# Multimodal fake news detection â€” complete project notebook
**Ali Abdulzahra | MSc project | Consolidated source and evidence companion**

This notebook brings together the project's data preparation, image audit and cleaning, unimodal training, fusion experiments, final holdout evaluation, explainability, later methodology checks and source-disjoint retraining. It includes the actual implementation rather than links to scripts alone.

The canonical code is the submission copy. Earlier local versions are retained in a labelled historical appendix. Consolidating the code does not mean the experiments were rerun: saved results are identified as saved evidence. The notebook was assembled with AI assistance from the existing project files; the report's AI-use section describes assistance during the project.

### How to use this notebook
1. **Read:** follow the sections in order; all Python source is visible.
2. **Run All for inspection:** cells beginning with `%%project_source` register source text without executing the experiment. The final checks compile that source and recompute the headline metrics from embedded saved predictions in a temporary folder. No GPU, original dataset or network is needed for these checks.
3. **Reproduce deliberately:** export a fresh working copy using the helper near the end, restore the external assets and choose individual scripts/stages. Training, downloads and analyses that write outputs are never automatically launched by Run All.

The inspection kernel needs Python, IPython and the standard library. Full experiments need their scientific/ML dependencies, data and weights. The embedded evidence supports inspection independently of the original F: drive; it does not include raw images or trained checkpoints.

### Contents
- [1. Research design and interpretation](#design)
- [2. Notebook machinery](#machinery)
- [3. Data preparation and cleaning](#data)
- [4. Unimodal baselines](#baselines)
- [5. Fusion experiments](#fusion)
- [6. Development diagnostics and explainability](#diagnostics)
- [7. Locked final holdout](#holdout)
- [8. Later methodology notebook](#methodology)
- [9. Source-disjoint retraining](#source)
- [10. Verification, configuration and historical sources](#support)
- [11. Saved evidence and reproduction controls](#reproduce)


<a id="design"></a>
## 1. Research design and interpretation

The research question is whether images add useful information to text for binary classification on cleaned Fakeddit samples. RoBERTa and ResNet-50 supply text and image baselines. Learned feature fusion and linear probes explore representations; probability fusion combines the two models' class-1 probabilities.

The image audit identified repeated regional-unavailability placeholders. Such files must be distinguished from valid duplicate content before filtering: a downloaded image can be readable yet semantically useless. Removal and failed-download patterns also affect which posts enter the multimodal subset. The code below records that selection rather than treating retained images as a random sample.

For late fusion, `p = alpha * p_text + (1 - alpha) * p_image`. Predictions are paired by post ID and checked for label agreement. Validation determines alpha; test data measures the frozen choice. Loading a test file before a search is different from using its labels in that search. The threshold is 0.50 for the ordinary locked evaluation.

The ordinary holdout has 5,000 cases and selects text weight 0.45 on development validation. Saved macro F1 is approximately 0.8000 (text), 0.7275 (image), and 0.8188 (fusion). The later source-disjoint experiment retrains on separate subreddit groups; its validation chooses text weight 0.00. On 2,739 test cases, macro F1 is approximately 0.7596 (text) and 0.6771 (image and locked fusion). Thus the ordinary gain does not establish reliable improvement on unseen sources.

The chronology is important: development results guided experiments; the ordinary frozen holdout is separate; later diagnostics and the source-disjoint experiment address further limitations. Creating a chronological manifest is not equivalent to training and evaluating a chronological model. Perceptual-hash matches are review candidates, not automatic proof of leakage. Fakeddit labels are dataset targets rather than independent fact-checking judgments.


<a id="machinery"></a>
## 2. Notebook machinery

The small cell magic below stores each source block under its original relative filename. Long files are split at top-level Python boundaries for readability and reassembled in order. Blank-line whitespace and line endings are normalised; Python statements are preserved. This preserves script entry points, command-line arguments, multiprocessing behaviour and separate namespaces. Editing a registered source block changes the exported working copy, not the original project. Restart and Run All after edits so the source registry is rebuilt consistently.

In [1]:
from pathlib import Path
import ast, base64, hashlib, io, json, os, subprocess, sys, tempfile, zipfile
from IPython.core.magic import register_cell_magic
from IPython.display import display, Markdown

SOURCE_PARTS = {}
@register_cell_magic
def project_source(line, cell):
    name, part = line.rsplit(" ", 1)
    SOURCE_PARTS.setdefault(name, {})[int(part)] = cell.rsplit("# END REGISTERED SOURCE BLOCK", 1)[0]

def registered_source(name):
    parts = SOURCE_PARTS[name]
    assert sorted(parts) == list(range(len(parts))), f"Missing source block: {name}"
    return "".join(parts[k] for k in sorted(parts))

print("Source registry ready. Experiment cells will be stored, not executed.")

Source registry ready. Experiment cells will be stored, not executed.


<a id="data"></a>
## 3. Data preparation and cleaning

Read the path constants and prerequisites before launching any stage. The ordering below follows the main dependencies; the code remains the authoritative record of each operation.

### 3.1 Audit fakeddit

Inspect dataset structure, labels, missing fields and sample counts before modelling.

**Source:** `multimodal-fake-news-detection/scripts/audit_fakeddit.py`  
**Imported modules:** `json`, `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/raw/fakeddit/multimodal_only_samples`
- `results/metrics`

The following cells contain the complete source; Run All registers it for inspection/export.

In [2]:
%%project_source multimodal-fake-news-detection/scripts/audit_fakeddit.py 0
from pathlib import Path
import json
import pandas as pd

BASE = Path("data/raw/fakeddit/multimodal_only_samples")

FILES = {
    "train": BASE / "multimodal_train.tsv",
    "validation": BASE / "multimodal_validate.tsv",
    "test": BASE / "multimodal_test_public.tsv",
}

OUTPUT_DIR = Path("results/metrics")
OUTPUT_DIR.mkdir(parents=True, exist_ok=True)

audit = {}

for split_name, path in FILES.items():
    print("=" * 80)
    print(f"{split_name.upper()}: {path}")
    print("=" * 80)

    df = pd.read_csv(path, sep="\t", low_memory=False)

    print(f"\nShape: {df.shape}")
    print(f"Memory: {df.memory_usage(deep=True).sum() / 1024**2:.2f} MB")

    print("\nColumns:")
    for column in df.columns:
        print(f"  - {column}")

    print("\nFirst 3 rows:")
    print(df.head(3).to_string())

    print("\nTop missing-value counts:")
    missing = df.isna().sum().sort_values(ascending=False)
    print(missing.head(20).to_string())

    print("\nLabel distributions:")
    label_info = {}

    for label_col in ["2_way_label", "3_way_label", "6_way_label"]:
        if label_col in df.columns:
            counts = df[label_col].value_counts(dropna=False).sort_index()
            print(f"\n{label_col}:")
            print(counts.to_string())

            label_info[label_col] = {
                str(k): int(v) for k, v in counts.items()
            }

    duplicate_info = {}

    for id_col in ["id", "submission_id"]:
        if id_col in df.columns:
            duplicate_info[id_col] = int(df[id_col].duplicated().sum())
            print(
                f"\nDuplicate {id_col} values: "
                f"{duplicate_info[id_col]}"
            )

    text_info = {}

    for text_col in ["clean_title", "title"]:
        if text_col in df.columns:
            lengths = df[text_col].fillna("").astype(str).str.len()

            text_info[text_col] = {
                "missing": int(df[text_col].isna().sum()),
                "empty": int((lengths == 0).sum()),
                "mean_length": float(lengths.mean()),
                "median_length": float(lengths.median()),
                "max_length": int(lengths.max()),
                "duplicates": int(df[text_col].duplicated().sum()),
            }

            print(f"\n{text_col} statistics:")
            for key, value in text_info[text_col].items():
                print(f"  {key}: {value}")

    image_info = {}

    for image_col in [
        "image_url",
        "hasImage",
        "image_id"
    ]:
        if image_col in df.columns:
            image_info[image_col] = {
                "missing": int(df[image_col].isna().sum()),
                "unique": int(df[image_col].nunique(dropna=True)),
            }

            print(f"\n{image_col}:")
            print(f"  missing: {image_info[image_col]['missing']}")
            print(f"  unique: {image_info[image_col]['unique']}")

    audit[split_name] = {
        "rows": int(len(df)),
        "columns": int(len(df.columns)),
        "column_names": list(df.columns),
        "memory_mb": float(
            df.memory_usage(deep=True).sum() / 1024**2
        ),
        "missing_values": {
            col: int(value)
            for col, value in missing.items()
        },
        "labels": label_info,
        "duplicates": duplicate_info,
        "text": text_info,
        "image": image_info,
    }

with open(
    OUTPUT_DIR / "fakeddit_audit.json",
    "w",
    encoding="utf-8"
) as f:
    json.dump(audit, f, indent=2)

print("\n" + "=" * 80)
print("Audit complete.")
print("Saved to results/metrics/fakeddit_audit.json")
print("=" * 80)
# END REGISTERED SOURCE BLOCK


### 3.2 Audit split leakage

Measure overlap across the official partitions before drawing independence conclusions.

**Source:** `multimodal-fake-news-detection/scripts/audit_split_leakage.py`  
**Imported modules:** `json`, `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/raw/fakeddit/multimodal_only_samples`
- `results/metrics/fakeddit_split_leakage.json`

The following cells contain the complete source; Run All registers it for inspection/export.

In [3]:
%%project_source multimodal-fake-news-detection/scripts/audit_split_leakage.py 0
from pathlib import Path
import json
import pandas as pd

BASE = Path("data/raw/fakeddit/multimodal_only_samples")

FILES = {
    "train": BASE / "multimodal_train.tsv",
    "validation": BASE / "multimodal_validate.tsv",
    "test": BASE / "multimodal_test_public.tsv",
}

OUTPUT = Path("results/metrics/fakeddit_split_leakage.json")
OUTPUT.parent.mkdir(parents=True, exist_ok=True)

USE_COLUMNS = [
    "id",
    "clean_title",
    "image_url",
    "2_way_label",
]

splits = {}

for name, path in FILES.items():
    print(f"Loading {name}...")
    splits[name] = pd.read_csv(
        path,
        sep="\t",
        usecols=USE_COLUMNS,
        low_memory=False
    )

pairs = [
    ("train", "validation"),
    ("train", "test"),
    ("validation", "test"),
]

report = {}

for left_name, right_name in pairs:
    left = splits[left_name]
    right = splits[right_name]

    print("\n" + "=" * 70)
    print(f"{left_name.upper()} vs {right_name.upper()}")
    print("=" * 70)

    pair_key = f"{left_name}_vs_{right_name}"
    report[pair_key] = {}

    # ID overlap
    left_ids = set(left["id"].dropna())
    right_ids = set(right["id"].dropna())
    id_overlap = left_ids.intersection(right_ids)

    print(f"ID overlap: {len(id_overlap)}")

    report[pair_key]["id_overlap"] = len(id_overlap)

    # Exact clean-title overlap
    left_titles = set(left["clean_title"].dropna())
    right_titles = set(right["clean_title"].dropna())
    title_overlap = left_titles.intersection(right_titles)

    print(f"Exact clean_title overlap: {len(title_overlap)}")

    report[pair_key]["clean_title_overlap"] = len(title_overlap)

    # Image URL overlap
    left_images = set(left["image_url"].dropna())
    right_images = set(right["image_url"].dropna())
    image_overlap = left_images.intersection(right_images)

    print(f"Image URL overlap: {len(image_overlap)}")

    report[pair_key]["image_url_overlap"] = len(image_overlap)

    # Exact text + image pair overlap
    left_pairs = set(
        zip(
            left["clean_title"].fillna(""),
            left["image_url"].fillna("")
        )
    )

    right_pairs = set(
        zip(
            right["clean_title"].fillna(""),
            right["image_url"].fillna("")
        )
    )

    pair_overlap = left_pairs.intersection(right_pairs)

    print(f"Exact text-image pair overlap: {len(pair_overlap)}")

    report[pair_key]["text_image_pair_overlap"] = len(pair_overlap)

with OUTPUT.open("w", encoding="utf-8") as f:
    json.dump(report, f, indent=2)

print("\nAudit complete.")
print(f"Saved to: {OUTPUT}")
# END REGISTERED SOURCE BLOCK


### 3.3 Prepare fakeddit

Read the release tables, standardise the fields and prepare processed splits, including the implemented duplicate-removal rules.

**Source:** `multimodal-fake-news-detection/scripts/prepare_fakeddit.py`  
**Imported modules:** `pandas`, `pathlib`  
**Top-level components:** `remove_training_duplicates`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/raw/fakeddit/multimodal_only_samples`
- `data/processed/fakeddit`

The following cells contain the complete source; Run All registers it for inspection/export.

In [4]:
%%project_source multimodal-fake-news-detection/scripts/prepare_fakeddit.py 0
from pathlib import Path
import pandas as pd

RAW = Path("data/raw/fakeddit/multimodal_only_samples")
OUT = Path("data/processed/fakeddit")
OUT.mkdir(parents=True, exist_ok=True)

FILES = {
    "train": RAW / "multimodal_train.tsv",
    "validation": RAW / "multimodal_validate.tsv",
    "test": RAW / "multimodal_test_public.tsv",
}

USECOLS = [
    "id",
    "clean_title",
    "image_url",
    "2_way_label",
]

processed = {}

for split, path in FILES.items():
    print(f"Processing {split}...")

    df = pd.read_csv(
        path,
        sep="\t",
        usecols=USECOLS,
        low_memory=False,
    )

    df = df.rename(
        columns={
            "clean_title": "text",
            "2_way_label": "label",
        }
    )

    df["split"] = split
    df["source_dataset"] = "fakeddit"

    df["text_length_chars"] = df["text"].str.len()
    df["text_length_words"] = (
        df["text"]
        .str.split()
        .str.len()
    )

    df["image_url_available"] = df["image_url"].notna()

    # Ensure expected types.
    df["id"] = df["id"].astype(str)
    df["text"] = df["text"].astype(str)
    df["label"] = df["label"].astype("int8")

    processed[split] = df

    print(f"  Rows: {len(df):,}")
    print(
        "  Labels:",
        df["label"].value_counts().sort_index().to_dict()
    )
    print(
        "  Missing image URLs:",
        int(df["image_url"].isna().sum())
    )

    df.to_parquet(
        OUT / f"{split}.parquet",
        index=False
    )

print("\nCreating leakage-reduced evaluation splits...")

train = processed["train"]
val = processed["validation"]
test = processed["test"]

train_titles = set(train["text"])
train_images = set(train["image_url"].dropna())

train_pairs = set(
    zip(
        train["text"],
        train["image_url"].fillna("")
    )
)

def remove_training_duplicates(df):
    pair_series = list(
        zip(
            df["text"],
            df["image_url"].fillna("")
        )
    )

    exact_pair_duplicate = pd.Series(
        [pair in train_pairs for pair in pair_series],
        index=df.index
    )

    cleaned = df.loc[~exact_pair_duplicate].copy()

    return cleaned, int(exact_pair_duplicate.sum())

val_clean, val_removed = remove_training_duplicates(val)
test_clean, test_removed = remove_training_duplicates(test)

val_clean.to_parquet(
    OUT / "validation_deduplicated.parquet",
    index=False
)

test_clean.to_parquet(
    OUT / "test_deduplicated.parquet",
    index=False
)

print(f"Validation exact pairs removed: {val_removed}")
print(f"Test exact pairs removed: {test_removed}")

print("\nProcessed files saved to:")
print(OUT)
# END REGISTERED SOURCE BLOCK


### 3.4 Create dev subset

Create the reproducible stratified development samples used for early experiments.

**Source:** `multimodal-fake-news-detection/scripts/create_dev_subset.py`  
**Imported modules:** `pandas`, `pathlib`, `sklearn`  
**Top-level components:** `stratified_sample`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit`
- `data/processed/fakeddit/development`

The following cells contain the complete source; Run All registers it for inspection/export.

In [5]:
%%project_source multimodal-fake-news-detection/scripts/create_dev_subset.py 0
from pathlib import Path

import pandas as pd
from sklearn.model_selection import train_test_split


SEED = 42

INPUT_DIR = Path("data/processed/fakeddit")
OUTPUT_DIR = Path("data/processed/fakeddit/development")

OUTPUT_DIR.mkdir(
    parents=True,
    exist_ok=True
)

TARGET_SIZES = {
    "train": 20_000,
    "validation": 3_000,
    "test": 3_000,
}

FILES = {
    "train": INPUT_DIR / "train.parquet",
    "validation": INPUT_DIR / "validation.parquet",
    "test": INPUT_DIR / "test.parquet",
}


def stratified_sample(df, sample_size):
    """
    Select a reproducible sample while preserving
    the binary label distribution.
    """

    if sample_size >= len(df):
        return df.copy()

    sampled, _ = train_test_split(
        df,
        train_size=sample_size,
        random_state=SEED,
        stratify=df["label"]
    )

    return (
        sampled
        .sample(frac=1, random_state=SEED)
        .reset_index(drop=True)
    )


for split_name, path in FILES.items():

    print("=" * 70)
    print(split_name.upper())
    print("=" * 70)

    df = pd.read_parquet(path)

    target_size = TARGET_SIZES[split_name]

    sampled = stratified_sample(
        df,
        target_size
    )

    original_distribution = (
        df["label"]
        .value_counts(normalize=True)
        .sort_index()
    )

    sampled_distribution = (
        sampled["label"]
        .value_counts(normalize=True)
        .sort_index()
    )

    print(f"Original size: {len(df):,}")
    print(f"Development size: {len(sampled):,}")

    print("\nOriginal label distribution:")
    print(original_distribution)

    print("\nDevelopment label distribution:")
    print(sampled_distribution)

    output_path = (
        OUTPUT_DIR /
        f"{split_name}.parquet"
    )

    sampled.to_parquet(
        output_path,
        index=False
    )

    print(f"\nSaved: {output_path}")

print("\nDevelopment subset complete.")
# END REGISTERED SOURCE BLOCK


### 3.5 Download dev images

Download development image candidates and record outcomes. This stage uses the network and writes images and logs.

**Source:** `multimodal-fake-news-detection/scripts/download_dev_images.py`  
**Imported modules:** `pandas`, `pathlib`, `requests`, `time`, `tqdm`  
**Top-level components:** `download_image`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development`
- `data/raw/fakeddit/development_images`
- `results/metrics`

The following cells contain the complete source; Run All registers it for inspection/export.

In [6]:
%%project_source multimodal-fake-news-detection/scripts/download_dev_images.py 0
from pathlib import Path
import time

import pandas as pd
import requests
from tqdm import tqdm


DATA_DIR = Path("data/processed/fakeddit/development")
IMAGE_ROOT = Path("data/raw/fakeddit/development_images")
LOG_DIR = Path("results/metrics")

IMAGE_ROOT.mkdir(parents=True, exist_ok=True)
LOG_DIR.mkdir(parents=True, exist_ok=True)

SPLITS = ["train", "validation", "test"]

TIMEOUT = 15
MAX_RETRIES = 3

HEADERS = {
    "User-Agent": (
        "Mozilla/5.0 "
        "(Windows NT 10.0; Win64; x64) "
        "AppleWebKit/537.36"
    )
}


def download_image(session, url, destination):
    """
    Download a single image with basic retry handling.
    """

    for attempt in range(1, MAX_RETRIES + 1):
        try:
            response = session.get(
                url,
                timeout=TIMEOUT,
                headers=HEADERS,
                stream=True
            )

            response.raise_for_status()

            content_type = response.headers.get(
                "Content-Type",
                ""
            ).lower()

            if "image" not in content_type:
                return False, f"non-image content: {content_type}"

            with destination.open("wb") as f:
                for chunk in response.iter_content(
                    chunk_size=8192
                ):
                    if chunk:
                        f.write(chunk)

            if destination.stat().st_size == 0:
                destination.unlink(missing_ok=True)
                return False, "zero-byte image"

            return True, ""

        except Exception as exc:
            if attempt == MAX_RETRIES:
                return False, str(exc)

            time.sleep(attempt * 1.5)

    return False, "unknown failure"


for split in SPLITS:

    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    manifest = pd.read_parquet(
        DATA_DIR / f"{split}.parquet"
    )

    image_dir = IMAGE_ROOT / split
    image_dir.mkdir(
        parents=True,
        exist_ok=True
    )

    failures = []
    skipped_missing_url = 0
    already_present = 0
    downloaded = 0

    with requests.Session() as session:

        for row in tqdm(
            manifest.itertuples(index=False),
            total=len(manifest),
            desc=f"Downloading {split}"
        ):

            sample_id = str(row.id)
            url = row.image_url

            destination = image_dir / f"{sample_id}.jpg"

            if destination.exists() and destination.stat().st_size > 0:
                already_present += 1
                continue

            if pd.isna(url) or not str(url).strip():
                skipped_missing_url += 1
                failures.append({
                    "id": sample_id,
                    "url": "",
                    "reason": "missing image URL"
                })
                continue

            success, reason = download_image(
                session,
                str(url),
                destination
            )

            if success:
                downloaded += 1
            else:
                destination.unlink(missing_ok=True)

                failures.append({
                    "id": sample_id,
                    "url": str(url),
                    "reason": reason
                })

    failure_df = pd.DataFrame(failures)

    failure_path = (
        LOG_DIR /
        f"fakeddit_{split}_image_download_failures.csv"
    )

    failure_df.to_csv(
        failure_path,
        index=False
    )

    print()
    print(f"Samples: {len(manifest):,}")
    print(f"Downloaded: {downloaded:,}")
    print(f"Already present: {already_present:,}")
    print(f"Missing URLs: {skipped_missing_url:,}")
    print(f"Failures: {len(failures):,}")
    print(f"Failure log: {failure_path}")

print("\nDevelopment image download complete.")
# END REGISTERED SOURCE BLOCK


### 3.6 Audit image integrity

Open downloaded images, calculate exact hashes and record unreadable or repeated files.

**Source:** `multimodal-fake-news-detection/scripts/audit_image_integrity.py`  
**Imported modules:** `PIL`, `hashlib`, `json`, `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/raw/fakeddit/development_images`
- `data/processed/fakeddit/development`
- `results/metrics`

The following cells contain the complete source; Run All registers it for inspection/export.

In [7]:
%%project_source multimodal-fake-news-detection/scripts/audit_image_integrity.py 0
from pathlib import Path
import hashlib
import json

import pandas as pd
from PIL import Image, UnidentifiedImageError


IMAGE_ROOT = Path("data/raw/fakeddit/development_images")
MANIFEST_ROOT = Path("data/processed/fakeddit/development")
OUTPUT_DIR = Path("results/metrics")
OUTPUT_DIR.mkdir(parents=True, exist_ok=True)

SPLITS = ["train", "validation", "test"]

summary = {}

for split in SPLITS:
    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    image_dir = IMAGE_ROOT / split
    manifest_path = MANIFEST_ROOT / f"{split}.parquet"

    manifest = pd.read_parquet(manifest_path)

    results = []
    hash_counts = {}

    for row in manifest.itertuples(index=False):
        sample_id = str(row.id)
        image_path = image_dir / f"{sample_id}.jpg"

        record = {
            "id": sample_id,
            "exists": image_path.exists(),
            "valid": False,
            "width": None,
            "height": None,
            "mode": None,
            "format": None,
            "size_bytes": None,
            "sha256": None,
            "error": None,
        }

        if not image_path.exists():
            record["error"] = "missing_file"
            results.append(record)
            continue

        try:
            record["size_bytes"] = image_path.stat().st_size

            with image_path.open("rb") as f:
                file_bytes = f.read()

            sha256 = hashlib.sha256(file_bytes).hexdigest()
            record["sha256"] = sha256

            hash_counts[sha256] = hash_counts.get(sha256, 0) + 1

            with Image.open(image_path) as img:
                img.verify()

            with Image.open(image_path) as img:
                img.load()

                record["width"] = img.width
                record["height"] = img.height
                record["mode"] = img.mode
                record["format"] = img.format

                if img.width <= 0 or img.height <= 0:
                    record["error"] = "invalid_dimensions"
                else:
                    record["valid"] = True

        except UnidentifiedImageError:
            record["error"] = "unidentified_image"

        except Exception as exc:
            record["error"] = str(exc)

        results.append(record)

    result_df = pd.DataFrame(results)

    duplicate_hashes = {
        h: count
        for h, count in hash_counts.items()
        if count > 1
    }

    output_csv = OUTPUT_DIR / f"fakeddit_{split}_image_integrity.csv"
    result_df.to_csv(output_csv, index=False)

    valid_count = int(result_df["valid"].sum())
    missing_count = int((~result_df["exists"]).sum())
    invalid_count = int(
        ((result_df["exists"]) & (~result_df["valid"])).sum()
    )

    suspicious_34641 = int(
        (result_df["size_bytes"] == 34641).sum()
    )

    duplicate_file_count = sum(
        count for count in duplicate_hashes.values()
    )

    print(f"Manifest rows: {len(result_df):,}")
    print(f"Valid images: {valid_count:,}")
    print(f"Missing files: {missing_count:,}")
    print(f"Invalid/corrupt images: {invalid_count:,}")
    print(f"Files exactly 34,641 bytes: {suspicious_34641:,}")
    print(f"Files involved in duplicate hashes: {duplicate_file_count:,}")
    print(f"Unique duplicated hashes: {len(duplicate_hashes):,}")

    summary[split] = {
        "manifest_rows": int(len(result_df)),
        "valid_images": valid_count,
        "missing_files": missing_count,
        "invalid_images": invalid_count,
        "files_34641_bytes": suspicious_34641,
        "duplicate_hash_groups": int(len(duplicate_hashes)),
        "files_in_duplicate_hash_groups": int(duplicate_file_count),
    }

with (OUTPUT_DIR / "fakeddit_image_integrity_summary.json").open(
    "w",
    encoding="utf-8"
) as f:
    json.dump(summary, f, indent=2)

print("\nImage integrity audit complete.")
# END REGISTERED SOURCE BLOCK


### 3.7 Inspect duplicate hashes

Inspect repeated image-hash groups to understand what the large duplicate group represents.

**Source:** `multimodal-fake-news-detection/scripts/inspect_duplicate_hashes.py`  
**Imported modules:** `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics`

The following cells contain the complete source; Run All registers it for inspection/export.

In [8]:
%%project_source multimodal-fake-news-detection/scripts/inspect_duplicate_hashes.py 0
from pathlib import Path
import pandas as pd

ROOT = Path("results/metrics")

for split in ["train", "validation", "test"]:
    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    path = ROOT / f"fakeddit_{split}_image_integrity.csv"
    df = pd.read_csv(path)

    valid = df[df["valid"] == True].copy()

    counts = (
        valid["sha256"]
        .value_counts()
        .reset_index()
    )

    counts.columns = ["sha256", "count"]

    repeated = counts[counts["count"] > 1]

    print("\nTop repeated hashes:")
    print(repeated.head(20).to_string(index=False))

    output = ROOT / f"fakeddit_{split}_duplicate_hashes.csv"
    repeated.to_csv(output, index=False)

    print(f"\nSaved: {output}")
# END REGISTERED SOURCE BLOCK


### 3.8 Create clean multimodal manifests

Build manifests for retained image/text pairs using the documented image-integrity exclusions.

**Source:** `multimodal-fake-news-detection/scripts/create_clean_multimodal_manifests.py`  
**Imported modules:** `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development`
- `results/metrics`
- `data/processed/fakeddit/development_clean`
- `data/raw/fakeddit/development_images`

The following cells contain the complete source; Run All registers it for inspection/export.

In [9]:
%%project_source multimodal-fake-news-detection/scripts/create_clean_multimodal_manifests.py 0
from pathlib import Path
import pandas as pd

MANIFEST_ROOT = Path("data/processed/fakeddit/development")
INTEGRITY_ROOT = Path("results/metrics")
OUTPUT_ROOT = Path("data/processed/fakeddit/development_clean")
OUTPUT_ROOT.mkdir(parents=True, exist_ok=True)

PLACEHOLDER_HASH = "faa24ec881e6040655c187a681d6dc496eb8aa41e1bd0652a180b3a40b457187"

for split in ["train", "validation", "test"]:
    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    manifest = pd.read_parquet(MANIFEST_ROOT / f"{split}.parquet")
    integrity = pd.read_csv(
        INTEGRITY_ROOT / f"fakeddit_{split}_image_integrity.csv"
    )

    integrity["id"] = integrity["id"].astype(str)
    manifest["id"] = manifest["id"].astype(str)

    integrity["is_placeholder"] = (
        integrity["sha256"] == PLACEHOLDER_HASH
    )

    integrity["image_usable"] = (
        integrity["exists"].eq(True)
        & integrity["valid"].eq(True)
        & ~integrity["is_placeholder"]
    )

    keep_cols = [
        "id",
        "exists",
        "valid",
        "image_usable",
        "is_placeholder",
        "width",
        "height",
        "size_bytes",
        "sha256",
        "error",
    ]

    merged = manifest.merge(
        integrity[keep_cols],
        on="id",
        how="left",
        validate="one_to_one"
    )

    merged["image_path"] = merged["id"].apply(
        lambda x: str(
            Path("data/raw/fakeddit/development_images")
            / split
            / f"{x}.jpg"
        )
    )

    usable = merged[merged["image_usable"] == True].copy()

    print(f"Original rows: {len(merged):,}")
    print(f"Usable multimodal rows: {len(usable):,}")
    print(f"Removed: {len(merged) - len(usable):,}")

    print("\nOriginal class distribution:")
    print(merged["label"].value_counts(normalize=True).sort_index())

    print("\nUsable class distribution:")
    print(usable["label"].value_counts(normalize=True).sort_index())

    merged.to_parquet(
        OUTPUT_ROOT / f"{split}_with_image_status.parquet",
        index=False
    )

    usable.to_parquet(
        OUTPUT_ROOT / f"{split}.parquet",
        index=False
    )

print("\nClean multimodal manifests complete.")
# END REGISTERED SOURCE BLOCK


### 3.9 Analyse placeholder sources

Examine the sources and labels associated with placeholder removals.

**Source:** `multimodal-fake-news-detection/scripts/analyse_placeholder_sources.py`  
**Imported modules:** `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/raw/fakeddit/multimodal_only_samples`
- `data/processed/fakeddit/development_clean`
- `results/metrics/fakeddit_placeholder_source_analysis.csv`

The following cells contain the complete source; Run All registers it for inspection/export.

In [10]:
%%project_source multimodal-fake-news-detection/scripts/analyse_placeholder_sources.py 0
from pathlib import Path
import pandas as pd

RAW_ROOT = Path("data/raw/fakeddit/multimodal_only_samples")
CLEAN_ROOT = Path("data/processed/fakeddit/development_clean")
OUTPUT = Path("results/metrics/fakeddit_placeholder_source_analysis.csv")

FILES = {
    "train": RAW_ROOT / "multimodal_train.tsv",
    "validation": RAW_ROOT / "multimodal_validate.tsv",
    "test": RAW_ROOT / "multimodal_test_public.tsv",
}

records = []

for split, raw_path in FILES.items():
    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    clean = pd.read_parquet(
        CLEAN_ROOT / f"{split}_with_image_status.parquet"
    )

    placeholder_ids = set(
        clean.loc[clean["is_placeholder"] == True, "id"].astype(str)
    )

    raw = pd.read_csv(
        raw_path,
        sep="\t",
        usecols=["id", "domain", "subreddit", "image_url"],
        low_memory=False
    )

    raw["id"] = raw["id"].astype(str)

    affected = raw[raw["id"].isin(placeholder_ids)].copy()

    print(f"Placeholder samples: {len(affected):,}")

    print("\nTop domains:")
    print(
        affected["domain"]
        .fillna("<missing>")
        .value_counts()
        .head(20)
        .to_string()
    )

    print("\nTop subreddits:")
    print(
        affected["subreddit"]
        .fillna("<missing>")
        .value_counts()
        .head(20)
        .to_string()
    )

    for domain, count in affected["domain"].fillna("<missing>").value_counts().items():
        records.append({
            "split": split,
            "domain": domain,
            "count": int(count)
        })

pd.DataFrame(records).to_csv(OUTPUT, index=False)

print(f"\nSaved: {OUTPUT}")
# END REGISTERED SOURCE BLOCK


### 3.10 Freeze fakeddit data

Record sample counts and ID fingerprints for the cleaned development partitions.

**Source:** `multimodal-fake-news-detection/scripts/freeze_fakeddit_data.py`  
**Imported modules:** `hashlib`, `json`, `pandas`, `pathlib`  
**Top-level components:** `hash_ids`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development_clean`
- `results/metrics/fakeddit_data_freeze.json`

The following cells contain the complete source; Run All registers it for inspection/export.

In [11]:
%%project_source multimodal-fake-news-detection/scripts/freeze_fakeddit_data.py 0
from pathlib import Path
import hashlib
import json

import pandas as pd


DATA_ROOT = Path("data/processed/fakeddit/development_clean")
OUTPUT = Path("results/metrics/fakeddit_data_freeze.json")

SPLITS = {
    "train": 13129,
    "validation": 1962,
    "test": 1965,
}


def hash_ids(ids):
    values = sorted(str(x) for x in ids)
    payload = "\n".join(values).encode("utf-8")
    return hashlib.sha256(payload).hexdigest()


summary = {}
id_sets = {}


for split, expected_count in SPLITS.items():

    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    path = DATA_ROOT / f"{split}.parquet"

    if not path.exists():
        raise FileNotFoundError(f"Missing dataset: {path}")

    df = pd.read_parquet(path)

    if len(df) != expected_count:
        raise ValueError(
            f"{split}: expected {expected_count:,} rows, "
            f"found {len(df):,}"
        )

    if df["id"].duplicated().any():
        raise ValueError(f"{split}: duplicate IDs detected.")

    labels = sorted(df["label"].unique().tolist())

    if labels != [0, 1]:
        raise ValueError(f"{split}: unexpected labels {labels}")

    if "image_usable" in df.columns:
        if not df["image_usable"].all():
            raise ValueError(f"{split}: unusable images remain.")

    missing_paths = 0

    if "image_path" in df.columns:
        missing_paths = sum(
            not Path(str(p)).exists()
            for p in df["image_path"]
        )

        if missing_paths:
            raise ValueError(
                f"{split}: {missing_paths} image paths do not exist."
            )

    ids = set(df["id"].astype(str))
    id_sets[split] = ids

    label_counts = (
        df["label"]
        .value_counts()
        .sort_index()
        .to_dict()
    )

    label_proportions = (
        df["label"]
        .value_counts(normalize=True)
        .sort_index()
        .to_dict()
    )

    split_hash = hash_ids(ids)

    summary[split] = {
        "rows": int(len(df)),
        "unique_ids": int(df["id"].nunique()),
        "label_counts": {
            str(k): int(v)
            for k, v in label_counts.items()
        },
        "label_proportions": {
            str(k): float(v)
            for k, v in label_proportions.items()
        },
        "sample_id_sha256": split_hash,
        "missing_image_paths": int(missing_paths),
    }

    print(f"Rows: {len(df):,}")
    print(f"Unique IDs: {df['id'].nunique():,}")
    print(f"Labels: {label_counts}")
    print(f"ID SHA256: {split_hash}")


train_val = id_sets["train"] & id_sets["validation"]
train_test = id_sets["train"] & id_sets["test"]
val_test = id_sets["validation"] & id_sets["test"]

summary["cross_split_id_overlap"] = {
    "train_validation": len(train_val),
    "train_test": len(train_test),
    "validation_test": len(val_test),
}

if train_val or train_test or val_test:
    raise ValueError("Cross-split ID overlap detected.")


OUTPUT.parent.mkdir(parents=True, exist_ok=True)

with OUTPUT.open("w", encoding="utf-8") as f:
    json.dump(summary, f, indent=2)

print("\n" + "=" * 70)
print("DATA FREEZE COMPLETE")
print("=" * 70)

print("\nCross-split ID overlap:")
print("Train / Validation:", len(train_val))
print("Train / Test:", len(train_test))
print("Validation / Test:", len(val_test))

print(f"\nFreeze record saved to: {OUTPUT}")
# END REGISTERED SOURCE BLOCK


### 3.11 Generate eda figures

Generate plots documenting dataset composition and image-cleaning effects.

**Source:** `multimodal-fake-news-detection/scripts/generate_eda_figures.py`  
**Imported modules:** `matplotlib`, `pandas`, `pathlib`  
**Top-level components:** `save_figure`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development`
- `data/processed/fakeddit/development_clean`
- `results/figures/eda`
- `results/metrics`

The following cells contain the complete source; Run All registers it for inspection/export.

In [12]:
%%project_source multimodal-fake-news-detection/scripts/generate_eda_figures.py 0
from pathlib import Path

import matplotlib.pyplot as plt
import pandas as pd


DEV_ROOT = Path("data/processed/fakeddit/development")
CLEAN_ROOT = Path("data/processed/fakeddit/development_clean")
FIGURE_ROOT = Path("results/figures/eda")
METRIC_ROOT = Path("results/metrics")

FIGURE_ROOT.mkdir(parents=True, exist_ok=True)
METRIC_ROOT.mkdir(parents=True, exist_ok=True)

SPLITS = ["train", "validation", "test"]

summary_rows = []


def save_figure(filename):
    plt.tight_layout()
    plt.savefig(FIGURE_ROOT / filename, dpi=300, bbox_inches="tight")
    plt.close()


# ============================================================
# Load datasets
# ============================================================

original = {}
status = {}
clean = {}

for split in SPLITS:
    original[split] = pd.read_parquet(
        DEV_ROOT / f"{split}.parquet"
    )

    status[split] = pd.read_parquet(
        CLEAN_ROOT / f"{split}_with_image_status.parquet"
    )

    clean[split] = pd.read_parquet(
        CLEAN_ROOT / f"{split}.parquet"
    )


# ============================================================
# 1. Original vs cleaned class distribution
# ============================================================

rows = []

for split in SPLITS:
    for dataset_name, df in [
        ("Original", original[split]),
        ("Cleaned", clean[split]),
    ]:
        counts = df["label"].value_counts().sort_index()

        for label, count in counts.items():
            rows.append({
                "split": split,
                "dataset": dataset_name,
                "label": int(label),
                "count": int(count),
                "proportion": count / len(df),
            })

class_df = pd.DataFrame(rows)

for split in SPLITS:
    subset = class_df[class_df["split"] == split]

    pivot = subset.pivot(
        index="label",
        columns="dataset",
        values="proportion"
    )

    ax = pivot.plot(kind="bar")

    ax.set_title(
        f"{split.capitalize()} class distribution: original vs cleaned"
    )
    ax.set_xlabel("Class label")
    ax.set_ylabel("Proportion")
    ax.set_ylim(0, 1)
    ax.legend(title="Dataset")

    plt.xticks(rotation=0)

    save_figure(
        f"{split}_class_distribution_original_vs_cleaned.png"
    )


# ============================================================
# 2. Image removal rate by class
# ============================================================

removal_rows = []

for split in SPLITS:
    df = status[split]

    removal = (
        df.groupby("label")["image_usable"]
        .apply(lambda x: 1 - x.mean())
    )

    for label, rate in removal.items():
        removal_rows.append({
            "split": split,
            "label": int(label),
            "removal_rate": float(rate),
        })

removal_df = pd.DataFrame(removal_rows)

pivot = removal_df.pivot(
    index="split",
    columns="label",
    values="removal_rate"
)

ax = pivot.plot(kind="bar")

ax.set_title("Unusable image rate by class and split")
ax.set_xlabel("Dataset split")
ax.set_ylabel("Removal rate")
ax.set_ylim(0, 1)
ax.legend(title="Class label")

plt.xticks(rotation=0)

save_figure("image_removal_rate_by_class.png")


# ============================================================
# 3. Overall usable image rate by split
# ============================================================

availability_rows = []

for split in SPLITS:
    df = status[split]

    usable = int(df["image_usable"].sum())
    total = len(df)

    availability_rows.append({
        "split": split,
        "usable": usable,
        "unusable": total - usable,
        "usable_rate": usable / total,
    })

availability_df = pd.DataFrame(availability_rows)

# END REGISTERED SOURCE BLOCK


In [13]:
%%project_source multimodal-fake-news-detection/scripts/generate_eda_figures.py 1
ax = availability_df.set_index("split")[
    ["usable", "unusable"]
].plot(
    kind="bar",
    stacked=True
)

ax.set_title("Usable and unusable images by split")
ax.set_xlabel("Dataset split")
ax.set_ylabel("Number of samples")

plt.xticks(rotation=0)

save_figure("usable_images_by_split.png")


# ============================================================
# 4. Text-length distribution
# ============================================================

combined_clean = pd.concat(
    [
        clean[split].assign(dataset_split=split)
        for split in SPLITS
    ],
    ignore_index=True
)

if "text_length_words" in combined_clean.columns:
    text_lengths = combined_clean["text_length_words"]
else:
    text_lengths = (
        combined_clean["text"]
        .fillna("")
        .astype(str)
        .str.split()
        .str.len()
    )

plt.figure()

plt.hist(
    text_lengths.clip(upper=text_lengths.quantile(0.995)),
    bins=50
)

plt.title("Text length distribution in cleaned multimodal dataset")
plt.xlabel("Number of words")
plt.ylabel("Number of samples")

save_figure("cleaned_text_length_distribution.png")


# ============================================================
# 5. Image width distribution
# ============================================================

image_rows = []

for split in SPLITS:
    df = status[split]

    usable = df[df["image_usable"] == True].copy()
    usable["dataset_split"] = split

    image_rows.append(usable)

usable_images = pd.concat(
    image_rows,
    ignore_index=True
)

width_limit = usable_images["width"].quantile(0.99)

plt.figure()

plt.hist(
    usable_images["width"].clip(upper=width_limit),
    bins=50
)

plt.title("Image width distribution")
plt.xlabel("Image width (pixels)")
plt.ylabel("Number of images")

save_figure("image_width_distribution.png")


# ============================================================
# 6. Image height distribution
# ============================================================

height_limit = usable_images["height"].quantile(0.99)

plt.figure()

plt.hist(
    usable_images["height"].clip(upper=height_limit),
    bins=50
)

plt.title("Image height distribution")
plt.xlabel("Image height (pixels)")
plt.ylabel("Number of images")

save_figure("image_height_distribution.png")


# ============================================================
# 7. Placeholder artefact counts
# ============================================================

placeholder_rows = []

for split in SPLITS:
    df = status[split]

    count = int(df["is_placeholder"].sum())

    placeholder_rows.append({
        "split": split,
        "placeholder_count": count,
    })

placeholder_df = pd.DataFrame(placeholder_rows)

ax = placeholder_df.set_index("split")[
    "placeholder_count"
].plot(kind="bar")

ax.set_title(
    "Repeated regional-unavailable placeholder images"
)
ax.set_xlabel("Dataset split")
ax.set_ylabel("Number of placeholder images")

plt.xticks(rotation=0)

save_figure("placeholder_images_by_split.png")


# ============================================================
# 8. Save numerical EDA summary
# ============================================================

for split in SPLITS:
    original_df = original[split]
    status_df = status[split]
    clean_df = clean[split]

    for label in sorted(original_df["label"].unique()):
        original_label = original_df[
            original_df["label"] == label
        ]

        status_label = status_df[
            status_df["label"] == label
        ]

        clean_label = clean_df[
            clean_df["label"] == label
        ]

        summary_rows.append({
            "split": split,
            "label": int(label),

            "original_count": len(original_label),
            "clean_count": len(clean_label),

            "original_proportion":
                len(original_label) / len(original_df),

            "clean_proportion":
                len(clean_label) / len(clean_df),

            "image_removal_rate":
                1 - status_label["image_usable"].mean(),

            "placeholder_count":
                int(status_label["is_placeholder"].sum()),
        })

# END REGISTERED SOURCE BLOCK


In [14]:
%%project_source multimodal-fake-news-detection/scripts/generate_eda_figures.py 2
summary_df = pd.DataFrame(summary_rows)

summary_df.to_csv(
    METRIC_ROOT / "fakeddit_eda_summary.csv",
    index=False
)


# ============================================================
# Console summary
# ============================================================

print("\n" + "=" * 70)
print("EDA COMPLETE")
print("=" * 70)

print("\nClean dataset sizes:")

for split in SPLITS:
    print(
        f"{split.capitalize():12s}: "
        f"{len(clean[split]):,}"
    )

print("\nFigures created:")

for figure in sorted(FIGURE_ROOT.glob("*.png")):
    print(f" - {figure}")

print(
    "\nSummary saved to:"
    "\nresults/metrics/fakeddit_eda_summary.csv"
)
# END REGISTERED SOURCE BLOCK


### 3.12 Audit token lengths

Measure token lengths to inform text truncation choices.

**Source:** `multimodal-fake-news-detection/scripts/audit_token_lengths.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `transformers`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit`
- `results/metrics/fakeddit_token_lengths.json`

The following cells contain the complete source; Run All registers it for inspection/export.

In [15]:
%%project_source multimodal-fake-news-detection/scripts/audit_token_lengths.py 0
from pathlib import Path
import json

import numpy as np
import pandas as pd
from transformers import AutoTokenizer


DATA_DIR = Path("data/processed/fakeddit")
OUTPUT = Path("results/metrics/fakeddit_token_lengths.json")

FILES = {
    "train": DATA_DIR / "train.parquet",
    "validation": DATA_DIR / "validation.parquet",
    "test": DATA_DIR / "test.parquet",
}

MODEL_NAME = "roberta-base"
BATCH_SIZE = 10000

print(f"Loading tokenizer: {MODEL_NAME}")

tokenizer = AutoTokenizer.from_pretrained(
    MODEL_NAME,
    use_fast=True
)

# Prevent warnings for long samples during the audit.
tokenizer.model_max_length = 1_000_000

report = {}

for split_name, path in FILES.items():

    print("\n" + "=" * 70)
    print(split_name.upper())
    print("=" * 70)

    df = pd.read_parquet(
        path,
        columns=["id", "text"]
    )

    lengths = []

    texts = df["text"].fillna("").astype(str).tolist()

    for start in range(0, len(texts), BATCH_SIZE):

        batch = texts[start:start + BATCH_SIZE]

        encoded = tokenizer(
            batch,
            add_special_tokens=True,
            padding=False,
            truncation=False,
            return_length=True
        )

        lengths.extend(encoded["length"])

        if start % 100000 == 0:
            print(
                f"Processed "
                f"{min(start + BATCH_SIZE, len(texts)):,}"
                f"/{len(texts):,}"
            )

    lengths = np.asarray(lengths)

    percentiles = {
        "p50": float(np.percentile(lengths, 50)),
        "p90": float(np.percentile(lengths, 90)),
        "p95": float(np.percentile(lengths, 95)),
        "p99": float(np.percentile(lengths, 99)),
        "p99_5": float(np.percentile(lengths, 99.5)),
        "p99_9": float(np.percentile(lengths, 99.9)),
    }

    thresholds = {}

    for threshold in [32, 64, 128, 256, 512]:
        percentage = (
            (lengths <= threshold).mean() * 100
        )

        thresholds[str(threshold)] = float(percentage)

    split_report = {
        "samples": int(len(lengths)),
        "mean": float(lengths.mean()),
        "median": float(np.median(lengths)),
        "min": int(lengths.min()),
        "max": int(lengths.max()),
        "percentiles": percentiles,
        "percentage_within_length": thresholds
    }

    report[split_name] = split_report

    print(f"Samples: {len(lengths):,}")
    print(f"Mean tokens: {lengths.mean():.2f}")
    print(f"Median tokens: {np.median(lengths):.0f}")
    print(f"Maximum tokens: {lengths.max()}")

    print("\nPercentiles:")

    for name, value in percentiles.items():
        print(f"  {name}: {value:.0f}")

    print("\nCoverage:")

    for threshold, percentage in thresholds.items():
        print(
            f"  <= {threshold:>3} tokens: "
            f"{percentage:.3f}%"
        )

OUTPUT.parent.mkdir(
    parents=True,
    exist_ok=True
)

with OUTPUT.open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        report,
        f,
        indent=2
    )

print("\n" + "=" * 70)
print("Token-length audit complete.")
print(f"Saved to: {OUTPUT}")
print("=" * 70)
# END REGISTERED SOURCE BLOCK


<a id="baselines"></a>
## 4. Unimodal baselines

Read the path constants and prerequisites before launching any stage. The ordering below follows the main dependencies; the code remains the authoritative record of each operation.

### 4.1 Train roberta baseline

Fine-tune the pretrained text encoder, evaluate validation performance and save the chosen checkpoint and metrics.

**Source:** `multimodal-fake-news-detection/scripts/train_roberta_baseline.py`  
**Imported modules:** `argparse`, `json`, `numpy`, `pandas`, `pathlib`, `random`, `sklearn`, `torch`, `transformers`  
**Top-level components:** `set_seed`, `TextDataset`, `compute_metrics`, `evaluate`, `train_epoch`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development_clean`
- `checkpoints/roberta_baseline`
- `results/metrics/roberta_baseline`

The following cells contain the complete source; Run All registers it for inspection/export.

In [16]:
%%project_source multimodal-fake-news-detection/scripts/train_roberta_baseline.py 0
import argparse
import json
import random
from pathlib import Path

import numpy as np
import pandas as pd
import torch

from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
    confusion_matrix,
)

from torch.optim import AdamW
from torch.utils.data import Dataset, DataLoader

from transformers import (
    AutoTokenizer,
    AutoModelForSequenceClassification,
    get_linear_schedule_with_warmup,
)


SEED = 42
MODEL_NAME = "roberta-base"
MAX_LENGTH = 64

DATA_ROOT = Path("data/processed/fakeddit/development_clean")
CHECKPOINT_ROOT = Path("checkpoints/roberta_baseline")
RESULT_ROOT = Path("results/metrics/roberta_baseline")

CHECKPOINT_ROOT.mkdir(parents=True, exist_ok=True)
RESULT_ROOT.mkdir(parents=True, exist_ok=True)


def set_seed(seed=SEED):
    random.seed(seed)
    np.random.seed(seed)

    torch.manual_seed(seed)

    if torch.cuda.is_available():
        torch.cuda.manual_seed_all(seed)

    torch.backends.cudnn.deterministic = True
    torch.backends.cudnn.benchmark = False


class TextDataset(Dataset):
    def __init__(self, dataframe, tokenizer):
        self.labels = torch.tensor(
            dataframe["label"].astype(int).values,
            dtype=torch.long
        )

        texts = (
            dataframe["text"]
            .fillna("")
            .astype(str)
            .tolist()
        )

        self.encodings = tokenizer(
            texts,
            padding="max_length",
            truncation=True,
            max_length=MAX_LENGTH,
            return_tensors="pt"
        )

    def __len__(self):
        return len(self.labels)

    def __getitem__(self, idx):
        item = {
            key: tensor[idx]
            for key, tensor in self.encodings.items()
        }

        item["labels"] = self.labels[idx]

        return item


def compute_metrics(labels, predictions, probabilities):
    metrics = {
        "accuracy": accuracy_score(labels, predictions),
        "precision": precision_score(
            labels,
            predictions,
            zero_division=0
        ),
        "recall": recall_score(
            labels,
            predictions,
            zero_division=0
        ),
        "f1": f1_score(
            labels,
            predictions,
            zero_division=0
        ),
        "f1_macro": f1_score(
        labels,
        predictions,
        average="macro",
        zero_division=0
        ),
    }

    try:
        metrics["roc_auc"] = roc_auc_score(
            labels,
            probabilities
        )
    except ValueError:
        metrics["roc_auc"] = None

    try:
        metrics["pr_auc"] = average_precision_score(
            labels,
            probabilities
        )
    except ValueError:
        metrics["pr_auc"] = None

    return metrics


def evaluate(model, loader, device):
    model.eval()

    total_loss = 0.0

    labels_all = []
    predictions_all = []
    probabilities_all = []

    with torch.no_grad():

        for batch in loader:

            labels = batch["labels"]

            batch = {
                key: value.to(device)
                for key, value in batch.items()
            }

            with torch.autocast(
                device_type="cuda",
                dtype=torch.float16,
                enabled=device.type == "cuda"
            ):
                outputs = model(**batch)

            loss = outputs.loss
            logits = outputs.logits

            total_loss += loss.item()

            probabilities = torch.softmax(
                logits,
                dim=1
            )[:, 1]

            predictions = torch.argmax(
                logits,
                dim=1
            )

            labels_all.extend(
                labels.cpu().numpy().tolist()
            )

            predictions_all.extend(
                predictions.cpu().numpy().tolist()
            )

            probabilities_all.extend(
                probabilities.cpu().numpy().tolist()
            )

    metrics = compute_metrics(
        labels_all,
        predictions_all,
        probabilities_all
    )

    metrics["loss"] = total_loss / len(loader)

    return (
        metrics,
        labels_all,
        predictions_all,
        probabilities_all
    )


# END REGISTERED SOURCE BLOCK


In [17]:
%%project_source multimodal-fake-news-detection/scripts/train_roberta_baseline.py 1
def train_epoch(
    model,
    loader,
    optimizer,
    scheduler,
    scaler,
    device
):
    model.train()

    total_loss = 0.0

    for step, batch in enumerate(loader, start=1):

        batch = {
            key: value.to(device)
            for key, value in batch.items()
        }

        optimizer.zero_grad(set_to_none=True)

        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=device.type == "cuda"
        ):
            outputs = model(**batch)
            loss = outputs.loss

        scaler.scale(loss).backward()

        scaler.unscale_(optimizer)

        torch.nn.utils.clip_grad_norm_(
            model.parameters(),
            max_norm=1.0
        )

        scaler.step(optimizer)
        scaler.update()

        scheduler.step()

        total_loss += loss.item()

        if step % 100 == 0:
            print(
                f"  Step {step:4d}/{len(loader)} "
                f"| Loss {total_loss / step:.4f}"
            )

    return total_loss / len(loader)


def main():

    parser = argparse.ArgumentParser()

    parser.add_argument(
        "--epochs",
        type=int,
        default=3
    )

    parser.add_argument(
        "--batch-size",
        type=int,
        default=16
    )

    parser.add_argument(
        "--lr",
        type=float,
        default=2e-5
    )

    parser.add_argument(
        "--smoke-test",
        action="store_true"
    )

    args = parser.parse_args()

    set_seed()

    device = torch.device(
        "cuda" if torch.cuda.is_available()
        else "cpu"
    )

    print("=" * 70)
    print("ROBERTA TEXT BASELINE")
    print("=" * 70)

    print(f"\nDevice: {device}")

    if device.type == "cuda":
        print(
            "GPU:",
            torch.cuda.get_device_name(0)
        )

    print(f"Model: {MODEL_NAME}")
    print(f"Max length: {MAX_LENGTH}")
    print(f"Batch size: {args.batch_size}")
    print(f"Learning rate: {args.lr}")
    print(f"Epochs: {args.epochs}")

    train_df = pd.read_parquet(
        DATA_ROOT / "train.parquet"
    )

    validation_df = pd.read_parquet(
        DATA_ROOT / "validation.parquet"
    )

    test_df = pd.read_parquet(
        DATA_ROOT / "test.parquet"
    )

    if args.smoke_test:

        print("\nSMOKE TEST MODE")

        train_df = train_df.sample(
            n=min(512, len(train_df)),
            random_state=SEED
        )

        validation_df = validation_df.sample(
            n=min(256, len(validation_df)),
            random_state=SEED
        )

        test_df = test_df.sample(
            n=min(256, len(test_df)),
            random_state=SEED
        )

        args.epochs = 1

    print("\nDataset sizes:")
    print(f"Train:      {len(train_df):,}")
    print(f"Validation: {len(validation_df):,}")
    print(f"Test:       {len(test_df):,}")

    tokenizer = AutoTokenizer.from_pretrained(
        MODEL_NAME
    )

    train_dataset = TextDataset(
        train_df,
        tokenizer
    )

    validation_dataset = TextDataset(
        validation_df,
        tokenizer
    )

    test_dataset = TextDataset(
        test_df,
        tokenizer
    )

    train_loader = DataLoader(
        train_dataset,
        batch_size=args.batch_size,
        shuffle=True,
        num_workers=0,
        pin_memory=device.type == "cuda"
    )

    validation_loader = DataLoader(
        validation_dataset,
        batch_size=args.batch_size,
        shuffle=False,
        num_workers=0,
        pin_memory=device.type == "cuda"
    )

    test_loader = DataLoader(
        test_dataset,
        batch_size=args.batch_size,
        shuffle=False,
        num_workers=0,
        pin_memory=device.type == "cuda"
    )

    model = AutoModelForSequenceClassification.from_pretrained(
        MODEL_NAME,
        num_labels=2
    )

    model.to(device)

    optimizer = AdamW(
        model.parameters(),
        lr=args.lr,
        weight_decay=0.01
    )

    total_steps = (
        len(train_loader)
        * args.epochs
    )

    warmup_steps = int(
        total_steps * 0.10
    )

    scheduler = get_linear_schedule_with_warmup(
        optimizer,
        num_warmup_steps=warmup_steps,
        num_training_steps=total_steps
    )

    scaler = torch.amp.GradScaler(
        "cuda",
        enabled=device.type == "cuda"
    )

    history = []

    best_f1 = -1.0
    epochs_without_improvement = 0
    patience = 2

    for epoch in range(
        1,
        args.epochs + 1
    ):

        print("\n" + "=" * 70)
        print(f"EPOCH {epoch}/{args.epochs}")
        print("=" * 70)

        train_loss = train_epoch(
            model,
            train_loader,
            optimizer,
            scheduler,
            scaler,
            device
        )

        val_metrics, _, _, _ = evaluate(
            model,
            validation_loader,
            device
        )

        print(
            f"\nTrain loss: {train_loss:.4f}"
        )

        print("\nValidation metrics:")

        for name, value in val_metrics.items():

            if value is None:
                print(f"{name:12s}: N/A")
            else:
                print(
                    f"{name:12s}: "
                    f"{value:.4f}"
                )

        epoch_record = {
            "epoch": epoch,
            "train_loss": train_loss,
            **{
                f"validation_{k}": v
                for k, v
                in val_metrics.items()
            }
        }

        history.append(epoch_record)

        current_f1 = val_metrics["f1_macro"]

        if current_f1 > best_f1:

            best_f1 = current_f1
            epochs_without_improvement = 0

            print(
                "\nNew best validation macro F1. "
                "Saving checkpoint."
            )

            model.save_pretrained(
                CHECKPOINT_ROOT
            )

            tokenizer.save_pretrained(
                CHECKPOINT_ROOT
            )

        else:

            epochs_without_improvement += 1

            print(
                "\nNo validation F1 improvement."
            )

            if (
                epochs_without_improvement
                >= patience
            ):

                print(
                    "Early stopping triggered."
                )

                break

    history_df = pd.DataFrame(history)

    history_df.to_csv(
        RESULT_ROOT / "training_history.csv",
        index=False
    )

    print("\nLoading best checkpoint...")

    best_model = (
        AutoModelForSequenceClassification
        .from_pretrained(
            CHECKPOINT_ROOT
        )
    )

    best_model.to(device)

    (
        test_metrics,
        test_labels,
        test_predictions,
        test_probabilities
    ) = evaluate(
        best_model,
        test_loader,
        device
    )

    print("\n" + "=" * 70)
    print("TEST RESULTS")
    print("=" * 70)

    for name, value in test_metrics.items():

        if value is None:
            print(f"{name:12s}: N/A")
        else:
            print(
                f"{name:12s}: "
                f"{value:.4f}"
            )

    matrix = confusion_matrix(
        test_labels,
        test_predictions
    )

    print("\nConfusion matrix:")
    print(matrix)

    with (
        RESULT_ROOT / "test_metrics.json"
    ).open(
        "w",
        encoding="utf-8"
    ) as f:

        json.dump(
            {
                **test_metrics,
                "confusion_matrix":
                    matrix.tolist(),
                "best_validation_f1":
                    best_f1,
                "model": MODEL_NAME,
                "max_length":
                    MAX_LENGTH,
                "seed":
                    SEED,
                "batch_size":
                    args.batch_size,
                "learning_rate":
                    args.lr,
            },
            f,
            indent=2
        )

    predictions_df = pd.DataFrame({
        "id": test_df["id"].astype(str),
        "label": test_labels,
        "prediction": test_predictions,
        "probability_class_1":
            test_probabilities
    })

    predictions_df.to_csv(
        RESULT_ROOT / "test_predictions.csv",
        index=False
    )

    print(
        "\nResults saved to:",
        RESULT_ROOT
    )

    print(
        "Best model saved to:",
        CHECKPOINT_ROOT
    )


# END REGISTERED SOURCE BLOCK


In [18]:
%%project_source multimodal-fake-news-detection/scripts/train_roberta_baseline.py 2
if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


### 4.2 Plot roberta baseline

Plot the stored text-model training/evaluation records.

**Source:** `multimodal-fake-news-detection/scripts/plot_roberta_baseline.py`  
**Imported modules:** `json`, `matplotlib`, `numpy`, `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/roberta_baseline`
- `results/figures/roberta_baseline`

The following cells contain the complete source; Run All registers it for inspection/export.

In [19]:
%%project_source multimodal-fake-news-detection/scripts/plot_roberta_baseline.py 0
from pathlib import Path

import json
import matplotlib.pyplot as plt
import pandas as pd
import numpy as np


RESULT_ROOT = Path("results/metrics/roberta_baseline")
FIGURE_ROOT = Path("results/figures/roberta_baseline")

FIGURE_ROOT.mkdir(parents=True, exist_ok=True)


# ------------------------------------------------------------
# Training history
# ------------------------------------------------------------

history = pd.read_csv(
    RESULT_ROOT / "training_history.csv"
)

plt.figure()

plt.plot(
    history["epoch"],
    history["train_loss"],
    marker="o",
    label="Training loss"
)

plt.plot(
    history["epoch"],
    history["validation_loss"],
    marker="o",
    label="Validation loss"
)

plt.xlabel("Epoch")
plt.ylabel("Loss")
plt.title("RoBERTa training and validation loss")
plt.xticks(history["epoch"])
plt.legend()

plt.tight_layout()
plt.savefig(
    FIGURE_ROOT / "training_validation_loss.png",
    dpi=300
)
plt.close()


# ------------------------------------------------------------
# Validation Macro F1
# ------------------------------------------------------------

plt.figure()

plt.plot(
    history["epoch"],
    history["validation_f1_macro"],
    marker="o"
)

plt.xlabel("Epoch")
plt.ylabel("Macro F1")
plt.title("RoBERTa validation Macro F1")
plt.xticks(history["epoch"])

plt.tight_layout()
plt.savefig(
    FIGURE_ROOT / "validation_macro_f1.png",
    dpi=300
)
plt.close()


# ------------------------------------------------------------
# Confusion matrix
# ------------------------------------------------------------

with (
    RESULT_ROOT / "test_metrics.json"
).open("r", encoding="utf-8") as f:
    metrics = json.load(f)

matrix = np.array(
    metrics["confusion_matrix"]
)

plt.figure()

plt.imshow(matrix)

plt.title("RoBERTa test confusion matrix")
plt.xlabel("Predicted class")
plt.ylabel("True class")

plt.xticks([0, 1], ["0", "1"])
plt.yticks([0, 1], ["0", "1"])

for i in range(2):
    for j in range(2):
        plt.text(
            j,
            i,
            str(matrix[i, j]),
            ha="center",
            va="center"
        )

plt.colorbar()

plt.tight_layout()
plt.savefig(
    FIGURE_ROOT / "test_confusion_matrix.png",
    dpi=300
)
plt.close()


print("RoBERTa baseline figures created.")

for path in sorted(FIGURE_ROOT.glob("*.png")):
    print(" -", path)
# END REGISTERED SOURCE BLOCK


### 4.3 Train resnet baseline

Train the image baseline on aligned clean samples and save checkpoints and evaluation records.

**Source:** `multimodal-fake-news-detection/scripts/train_resnet_baseline.py`  
**Imported modules:** `PIL`, `argparse`, `json`, `numpy`, `pandas`, `pathlib`, `random`, `sklearn`, `torch`, `torchvision`  
**Top-level components:** `set_seed`, `ImageDataset`, `compute_metrics`, `evaluate`, `train_epoch`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development_clean`
- `checkpoints/resnet50_baseline`
- `results/metrics/resnet50_baseline`

The following cells contain the complete source; Run All registers it for inspection/export.

In [20]:
%%project_source multimodal-fake-news-detection/scripts/train_resnet_baseline.py 0
import argparse
import json
import random
from pathlib import Path

import numpy as np
import pandas as pd
from PIL import Image

import torch
import torch.nn as nn

from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
    confusion_matrix,
)

from torch.optim import AdamW
from torch.utils.data import Dataset, DataLoader

from torchvision.models import (
    resnet50,
    ResNet50_Weights,
)

from torchvision import transforms


SEED = 42

DATA_ROOT = Path("data/processed/fakeddit/development_clean")
CHECKPOINT_ROOT = Path("checkpoints/resnet50_baseline")
RESULT_ROOT = Path("results/metrics/resnet50_baseline")

CHECKPOINT_ROOT.mkdir(parents=True, exist_ok=True)
RESULT_ROOT.mkdir(parents=True, exist_ok=True)


def set_seed(seed=SEED):
    random.seed(seed)
    np.random.seed(seed)

    torch.manual_seed(seed)

    if torch.cuda.is_available():
        torch.cuda.manual_seed_all(seed)

    torch.backends.cudnn.deterministic = True
    torch.backends.cudnn.benchmark = False


class ImageDataset(Dataset):
    def __init__(self, dataframe, transform):
        self.df = dataframe.reset_index(drop=True)
        self.transform = transform

    def __len__(self):
        return len(self.df)

    def __getitem__(self, idx):

        row = self.df.iloc[idx]

        image_path = Path(str(row["image_path"]))

        with Image.open(image_path) as image:
            image = image.convert("RGB")

        image = self.transform(image)

        label = torch.tensor(
            int(row["label"]),
            dtype=torch.long
        )

        return {
            "image": image,
            "label": label
        }


def compute_metrics(
    labels,
    predictions,
    probabilities
):
    metrics = {
        "accuracy": accuracy_score(
            labels,
            predictions
        ),

        "precision": precision_score(
            labels,
            predictions,
            zero_division=0
        ),

        "recall": recall_score(
            labels,
            predictions,
            zero_division=0
        ),

        "f1": f1_score(
            labels,
            predictions,
            zero_division=0
        ),

        "f1_macro": f1_score(
            labels,
            predictions,
            average="macro",
            zero_division=0
        ),
    }

    try:
        metrics["roc_auc"] = roc_auc_score(
            labels,
            probabilities
        )
    except ValueError:
        metrics["roc_auc"] = None

    try:
        metrics["pr_auc"] = average_precision_score(
            labels,
            probabilities
        )
    except ValueError:
        metrics["pr_auc"] = None

    return metrics


def evaluate(
    model,
    loader,
    device
):
    model.eval()

    total_loss = 0.0

    labels_all = []
    predictions_all = []
    probabilities_all = []

    criterion = nn.CrossEntropyLoss()

    with torch.no_grad():

        for batch in loader:

            images = batch["image"].to(
                device,
                non_blocking=True
            )

            labels = batch["label"].to(
                device,
                non_blocking=True
            )

            with torch.autocast(
                device_type="cuda",
                dtype=torch.float16,
                enabled=device.type == "cuda"
            ):

                logits = model(images)

                loss = criterion(
                    logits,
                    labels
                )

            probabilities = torch.softmax(
                logits,
                dim=1
            )[:, 1]

            predictions = torch.argmax(
                logits,
                dim=1
            )

            total_loss += loss.item()

            labels_all.extend(
                labels.cpu().numpy().tolist()
            )

            predictions_all.extend(
                predictions.cpu().numpy().tolist()
            )

            probabilities_all.extend(
                probabilities.cpu().numpy().tolist()
            )

    metrics = compute_metrics(
        labels_all,
        predictions_all,
        probabilities_all
    )

    metrics["loss"] = (
        total_loss / len(loader)
    )

    return (
        metrics,
        labels_all,
        predictions_all,
        probabilities_all
    )


# END REGISTERED SOURCE BLOCK


In [21]:
%%project_source multimodal-fake-news-detection/scripts/train_resnet_baseline.py 1
def train_epoch(
    model,
    loader,
    optimizer,
    scaler,
    criterion,
    device
):
    model.train()

    total_loss = 0.0

    for step, batch in enumerate(
        loader,
        start=1
    ):

        images = batch["image"].to(
            device,
            non_blocking=True
        )

        labels = batch["label"].to(
            device,
            non_blocking=True
        )

        optimizer.zero_grad(
            set_to_none=True
        )

        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=device.type == "cuda"
        ):

            logits = model(images)

            loss = criterion(
                logits,
                labels
            )

        scaler.scale(loss).backward()

        scaler.unscale_(
            optimizer
        )

        torch.nn.utils.clip_grad_norm_(
            model.parameters(),
            max_norm=1.0
        )

        scaler.step(
            optimizer
        )

        scaler.update()

        total_loss += loss.item()

        if step % 100 == 0:

            print(
                f"  Step {step:4d}/{len(loader)} "
                f"| Loss {total_loss / step:.4f}"
            )

    return (
        total_loss / len(loader)
    )


def main():

    parser = argparse.ArgumentParser()

    parser.add_argument(
        "--epochs",
        type=int,
        default=3
    )

    parser.add_argument(
        "--batch-size",
        type=int,
        default=32
    )

    parser.add_argument(
        "--lr",
        type=float,
        default=1e-4
    )

    parser.add_argument(
        "--num-workers",
        type=int,
        default=4
    )

    parser.add_argument(
        "--smoke-test",
        action="store_true"
    )

    args = parser.parse_args()

    set_seed()

    device = torch.device(
        "cuda"
        if torch.cuda.is_available()
        else "cpu"
    )

    if args.smoke_test:
        args.epochs = 1

    print("=" * 70)
    print("RESNET-50 IMAGE BASELINE")
    print("=" * 70)

    print(f"\nDevice: {device}")

    if device.type == "cuda":
        print(
            "GPU:",
            torch.cuda.get_device_name(0)
        )

    print("Model: ResNet-50")
    print("Input size: 224 x 224")
    print(f"Batch size: {args.batch_size}")
    print(f"Learning rate: {args.lr}")
    print(f"Epochs: {args.epochs}")
    print(
        f"DataLoader workers: "
        f"{args.num_workers}"
    )

    train_df = pd.read_parquet(
        DATA_ROOT / "train.parquet"
    )

    validation_df = pd.read_parquet(
        DATA_ROOT / "validation.parquet"
    )

    test_df = pd.read_parquet(
        DATA_ROOT / "test.parquet"
    )

    if args.smoke_test:

        print("\nSMOKE TEST MODE")

        train_df = train_df.sample(
            n=min(512, len(train_df)),
            random_state=SEED
        )

        validation_df = validation_df.sample(
            n=min(256, len(validation_df)),
            random_state=SEED
        )

        test_df = test_df.sample(
            n=min(256, len(test_df)),
            random_state=SEED
        )

    print("\nDataset sizes:")

    print(
        f"Train:      {len(train_df):,}"
    )

    print(
        f"Validation: {len(validation_df):,}"
    )

    print(
        f"Test:       {len(test_df):,}"
    )


    # --------------------------------------------------------
    # Image preprocessing
    # --------------------------------------------------------

    transform = transforms.Compose([
        transforms.Resize(
            (224, 224)
        ),

        transforms.ToTensor(),

        transforms.Normalize(
            mean=[
                0.485,
                0.456,
                0.406
            ],
            std=[
                0.229,
                0.224,
                0.225
            ]
        ),
    ])


    train_dataset = ImageDataset(
        train_df,
        transform
    )

    validation_dataset = ImageDataset(
        validation_df,
        transform
    )

    test_dataset = ImageDataset(
        test_df,
        transform
    )


    loader_kwargs = {
        "num_workers":
            args.num_workers,

        "pin_memory":
            device.type == "cuda",
    }

    if args.num_workers > 0:
        loader_kwargs[
            "persistent_workers"
        ] = True


    train_loader = DataLoader(
        train_dataset,
        batch_size=args.batch_size,
        shuffle=True,
        **loader_kwargs
    )

    validation_loader = DataLoader(
        validation_dataset,
        batch_size=args.batch_size,
        shuffle=False,
        **loader_kwargs
    )

    test_loader = DataLoader(
        test_dataset,
        batch_size=args.batch_size,
        shuffle=False,
        **loader_kwargs
    )


    # --------------------------------------------------------
    # Pretrained ResNet
    # --------------------------------------------------------

    weights = (
        ResNet50_Weights.IMAGENET1K_V2
    )

    model = resnet50(
        weights=weights
    )

    num_features = (
        model.fc.in_features
    )

    model.fc = nn.Linear(
        num_features,
        2
    )

    model.to(device)


    criterion = (
        nn.CrossEntropyLoss()
    )


    optimizer = AdamW(
        model.parameters(),
        lr=args.lr,
        weight_decay=0.01
    )


    scaler = torch.amp.GradScaler(
        "cuda",
        enabled=device.type == "cuda"
    )


    history = []

    best_macro_f1 = -1.0
    epochs_without_improvement = 0

    patience = 2


    # --------------------------------------------------------
    # Training
    # --------------------------------------------------------

    for epoch in range(
        1,
        args.epochs + 1
    ):

        print("\n" + "=" * 70)

        print(
            f"EPOCH {epoch}/{args.epochs}"
        )

        print("=" * 70)


        train_loss = train_epoch(
            model,
            train_loader,
            optimizer,
            scaler,
            criterion,
            device
        )


        (
            val_metrics,
            _,
            _,
            _
        ) = evaluate(
            model,
            validation_loader,
            device
        )


        print(
            f"\nTrain loss: "
            f"{train_loss:.4f}"
        )


        print(
            "\nValidation metrics:"
        )


        for name, value in (
            val_metrics.items()
        ):

            if value is None:

                print(
                    f"{name:12s}: N/A"
                )

            else:

                print(
                    f"{name:12s}: "
                    f"{value:.4f}"
                )


        history.append({
            "epoch": epoch,
            "train_loss": train_loss,

            **{
                f"validation_{key}":
                    value

                for key, value
                in val_metrics.items()
            }
        })


        current_macro_f1 = (
            val_metrics["f1_macro"]
        )


        if (
            current_macro_f1
            > best_macro_f1
        ):

            best_macro_f1 = (
                current_macro_f1
            )

            epochs_without_improvement = 0


            print(
                "\nNew best validation "
                "macro F1. "
                "Saving checkpoint."
            )


            torch.save(
                {
                    "model_state_dict":
                        model.state_dict(),

                    "model":
                        "resnet50",

                    "num_classes":
                        2,

                    "validation_macro_f1":
                        best_macro_f1,
                },

                CHECKPOINT_ROOT
                / "best_model.pt"
            )


        else:

            epochs_without_improvement += 1

            print(
                "\nNo validation macro "
                "F1 improvement."
            )


            if (
                epochs_without_improvement
                >= patience
            ):

                print(
                    "Early stopping "
                    "triggered."
                )

                break


    # --------------------------------------------------------
    # Save training history
    # --------------------------------------------------------

    pd.DataFrame(
        history
    ).to_csv(
        RESULT_ROOT
        / "training_history.csv",
        index=False
    )


    # --------------------------------------------------------
    # Load best checkpoint
    # --------------------------------------------------------

    print(
        "\nLoading best checkpoint..."
    )


    checkpoint = torch.load(
        CHECKPOINT_ROOT
        / "best_model.pt",
        map_location=device,
        weights_only=True
    )


    model.load_state_dict(
        checkpoint[
            "model_state_dict"
        ]
    )


    # --------------------------------------------------------
    # Final test evaluation
    # --------------------------------------------------------

    (
        test_metrics,
        test_labels,
        test_predictions,
        test_probabilities
    ) = evaluate(
        model,
        test_loader,
        device
    )


    print("\n" + "=" * 70)
    print("TEST RESULTS")
    print("=" * 70)


    for name, value in (
        test_metrics.items()
    ):

        if value is None:

            print(
                f"{name:12s}: N/A"
            )

        else:

            print(
                f"{name:12s}: "
                f"{value:.4f}"
            )


    matrix = confusion_matrix(
        test_labels,
        test_predictions
    )


    print(
        "\nConfusion matrix:"
    )

    print(matrix)


    # --------------------------------------------------------
    # Save metrics
    # --------------------------------------------------------

    with (
        RESULT_ROOT
        / "test_metrics.json"
    ).open(
        "w",
        encoding="utf-8"
    ) as f:

        json.dump(
            {
                **test_metrics,

                "confusion_matrix":
                    matrix.tolist(),

                "best_validation_macro_f1":
                    best_macro_f1,

                "model":
                    "resnet50",

                "weights":
                    "IMAGENET1K_V2",

                "image_size":
                    224,

                "seed":
                    SEED,

                "batch_size":
                    args.batch_size,

                "learning_rate":
                    args.lr,
            },

            f,
            indent=2
        )


    predictions_df = pd.DataFrame({
        "id":
            test_df["id"].astype(str),

        "label":
            test_labels,

        "prediction":
            test_predictions,

        "probability_class_1":
            test_probabilities
    })


    predictions_df.to_csv(
        RESULT_ROOT
        / "test_predictions.csv",
        index=False
    )


    print(
        "\nResults saved to:",
        RESULT_ROOT
    )

    print(
        "Best model saved to:",
        CHECKPOINT_ROOT
    )


# END REGISTERED SOURCE BLOCK


In [22]:
%%project_source multimodal-fake-news-detection/scripts/train_resnet_baseline.py 2
if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


<a id="fusion"></a>
## 5. Fusion experiments

Feature fusion consumes exported representations; probability fusion consumes per-ID probabilities. Training or tuning a fusion head is not interchangeable with selecting the late-fusion coefficient.

### 5.1 Extract multimodal features

Use trained encoders to export aligned text and image representations for fusion experiments.

**Source:** `multimodal-fake-news-detection/scripts/extract_multimodal_features.py`  
**Imported modules:** `PIL`, `argparse`, `pandas`, `pathlib`, `torch`, `torchvision`, `transformers`  
**Top-level components:** `MultimodalDataset`, `load_roberta`, `load_resnet`, `extract_split`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development_clean`
- `checkpoints/roberta_baseline`
- `checkpoints/resnet50_baseline/best_model.pt`
- `data/processed/fakeddit/multimodal_features`
- `data/processed/fakeddit/multimodal_features_smoke`

The following cells contain the complete source; Run All registers it for inspection/export.

In [23]:
%%project_source multimodal-fake-news-detection/scripts/extract_multimodal_features.py 0
import argparse
from pathlib import Path

import pandas as pd
from PIL import Image

import torch
import torch.nn as nn
from torch.utils.data import Dataset, DataLoader

from transformers import (
    AutoTokenizer,
    AutoModelForSequenceClassification,
)

from torchvision.models import resnet50
from torchvision import transforms


SEED = 42
MAX_LENGTH = 64

DATA_ROOT = Path("data/processed/fakeddit/development_clean")

ROBERTA_CHECKPOINT = Path("checkpoints/roberta_baseline")
RESNET_CHECKPOINT = Path("checkpoints/resnet50_baseline/best_model.pt")

OUTPUT_ROOT = Path("data/processed/fakeddit/multimodal_features")


class MultimodalDataset(Dataset):

    def __init__(
        self,
        dataframe,
        tokenizer,
        image_transform
    ):
        self.df = dataframe.reset_index(drop=True)

        self.tokenizer = tokenizer
        self.image_transform = image_transform

    def __len__(self):
        return len(self.df)

    def __getitem__(self, idx):

        row = self.df.iloc[idx]

        sample_id = str(row["id"])

        text = str(row["text"])

        tokens = self.tokenizer(
            text,
            truncation=True,
            max_length=MAX_LENGTH,
            padding="max_length",
            return_tensors="pt"
        )

        tokens = {
            key: value.squeeze(0)
            for key, value in tokens.items()
        }

        image_path = Path(
            str(row["image_path"])
        )

        with Image.open(image_path) as image:
            image = image.convert("RGB")
            image = self.image_transform(image)

        label = int(row["label"])

        return {
            "id": sample_id,
            "input_ids": tokens["input_ids"],
            "attention_mask": tokens["attention_mask"],
            "image": image,
            "label": label,
        }


def load_roberta(device):

    print("Loading fine-tuned RoBERTa...")

    model = (
        AutoModelForSequenceClassification
        .from_pretrained(
            ROBERTA_CHECKPOINT
        )
    )

    model.to(device)
    model.eval()

    for parameter in model.parameters():
        parameter.requires_grad = False

    return model


def load_resnet(device):

    print("Loading fine-tuned ResNet-50...")

    checkpoint = torch.load(
        RESNET_CHECKPOINT,
        map_location="cpu",
        weights_only=True
    )

    model = resnet50(
        weights=None
    )

    num_features = model.fc.in_features

    model.fc = nn.Linear(
        num_features,
        2
    )

    model.load_state_dict(
        checkpoint["model_state_dict"]
    )

    # Remove classifier so output becomes
    # the 2048-dimensional visual feature vector.
    model.fc = nn.Identity()

    model.to(device)
    model.eval()

    for parameter in model.parameters():
        parameter.requires_grad = False

    return model


@torch.no_grad()
def extract_split(
    split,
    dataframe,
    tokenizer,
    roberta,
    resnet,
    image_transform,
    device,
    batch_size,
    num_workers,
    output_root
):

    print("\n" + "=" * 70)
    print(split.upper())
    print("=" * 70)

    dataset = MultimodalDataset(
        dataframe,
        tokenizer,
        image_transform
    )

    loader_kwargs = {
        "batch_size": batch_size,
        "shuffle": False,
        "num_workers": num_workers,
        "pin_memory": device.type == "cuda",
    }

    if num_workers > 0:
        loader_kwargs[
            "persistent_workers"
        ] = True

    loader = DataLoader(
        dataset,
        **loader_kwargs
    )

    all_ids = []
    all_labels = []

    all_text_features = []
    all_image_features = []

    for step, batch in enumerate(
        loader,
        start=1
    ):

        input_ids = batch[
            "input_ids"
        ].to(
            device,
            non_blocking=True
        )

        attention_mask = batch[
            "attention_mask"
        ].to(
            device,
            non_blocking=True
        )

        images = batch[
            "image"
        ].to(
            device,
            non_blocking=True
        )

        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=device.type == "cuda"
        ):

            roberta_output = (
                roberta.roberta(
                    input_ids=input_ids,
                    attention_mask=attention_mask
                )
            )

            # First-token representation
            text_features = (
                roberta_output
                .last_hidden_state[:, 0, :]
            )

            image_features = resnet(
                images
            )

        all_text_features.append(
            text_features.float().cpu()
        )

        all_image_features.append(
            image_features.float().cpu()
        )

        all_labels.append(
            batch["label"].long()
        )

        all_ids.extend(
            batch["id"]
        )

        if step % 100 == 0:
            print(
                f"  Batch {step:4d}/{len(loader)}"
            )

    text_features = torch.cat(
        all_text_features,
        dim=0
    )

    image_features = torch.cat(
        all_image_features,
        dim=0
    )

    labels = torch.cat(
        all_labels,
        dim=0
    )

    if text_features.shape[0] != len(dataframe):
        raise ValueError(
            "Text feature row count mismatch."
        )

    if image_features.shape[0] != len(dataframe):
        raise ValueError(
            "Image feature row count mismatch."
        )

    print(
        f"\nSamples:        {len(all_ids):,}"
    )

    print(
        "Text features: ",
        tuple(text_features.shape)
    )

    print(
        "Image features:",
        tuple(image_features.shape)
    )

    output_root.mkdir(
        parents=True,
        exist_ok=True
    )

    output_path = (
        output_root
        / f"{split}.pt"
    )

    torch.save(
        {
            "ids": all_ids,
            "labels": labels,
            "text_features":
                text_features,
            "image_features":
                image_features,
        },
        output_path
    )

    print(
        f"Saved: {output_path}"
    )


# END REGISTERED SOURCE BLOCK


In [24]:
%%project_source multimodal-fake-news-detection/scripts/extract_multimodal_features.py 1
def main():

    parser = argparse.ArgumentParser()

    parser.add_argument(
        "--batch-size",
        type=int,
        default=32
    )

    parser.add_argument(
        "--num-workers",
        type=int,
        default=4
    )

    parser.add_argument(
        "--smoke-test",
        action="store_true"
    )

    args = parser.parse_args()

    torch.manual_seed(SEED)

    device = torch.device(
        "cuda"
        if torch.cuda.is_available()
        else "cpu"
    )

    print("=" * 70)
    print("MULTIMODAL FEATURE EXTRACTION")
    print("=" * 70)

    print(f"\nDevice: {device}")

    if device.type == "cuda":
        print(
            "GPU:",
            torch.cuda.get_device_name(0)
        )

    tokenizer = (
        AutoTokenizer
        .from_pretrained(
            ROBERTA_CHECKPOINT
        )
    )

    roberta = load_roberta(
        device
    )

    resnet = load_resnet(
        device
    )

    image_transform = transforms.Compose([
        transforms.Resize(
            (224, 224)
        ),

        transforms.ToTensor(),

        transforms.Normalize(
            mean=[
                0.485,
                0.456,
                0.406
            ],
            std=[
                0.229,
                0.224,
                0.225
            ]
        ),
    ])

    output_root = OUTPUT_ROOT

    if args.smoke_test:

        print("\nSMOKE TEST MODE")

        output_root = Path(
            "data/processed/fakeddit/"
            "multimodal_features_smoke"
        )

    for split in [
        "train",
        "validation",
        "test"
    ]:

        df = pd.read_parquet(
            DATA_ROOT / f"{split}.parquet"
        )

        if args.smoke_test:

            df = df.sample(
                n=min(256, len(df)),
                random_state=SEED
            ).reset_index(drop=True)

        extract_split(
            split=split,
            dataframe=df,
            tokenizer=tokenizer,
            roberta=roberta,
            resnet=resnet,
            image_transform=image_transform,
            device=device,
            batch_size=args.batch_size,
            num_workers=args.num_workers,
            output_root=output_root
        )

    print("\n" + "=" * 70)
    print("FEATURE EXTRACTION COMPLETE")
    print("=" * 70)


if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


### 5.2 Train multimodal fusion

Train a fusion MLP on extracted representations, including the implemented standardisation and regularisation controls.

**Source:** `multimodal-fake-news-detection/scripts/train_multimodal_fusion.py`  
**Imported modules:** `argparse`, `json`, `numpy`, `pandas`, `pathlib`, `random`, `sklearn`, `torch`  
**Top-level components:** `set_seed`, `load_features`, `standardize`, `FusionMLP`, `compute_metrics`, `evaluate`, `train_epoch`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/multimodal_features`
- `checkpoints/multimodal_fusion_baseline`
- `results/metrics/multimodal_fusion_baseline`

The following cells contain the complete source; Run All registers it for inspection/export.

In [25]:
%%project_source multimodal-fake-news-detection/scripts/train_multimodal_fusion.py 0
import argparse
import json
import random
from pathlib import Path

import numpy as np
import pandas as pd
import torch
import torch.nn as nn

from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
    confusion_matrix,
)

from torch.optim import AdamW
from torch.utils.data import TensorDataset, DataLoader


SEED = 42

FEATURE_ROOT = Path(
    "data/processed/fakeddit/multimodal_features"
)

CHECKPOINT_ROOT = Path(
    "checkpoints/multimodal_fusion_baseline"
)

RESULT_ROOT = Path(
    "results/metrics/multimodal_fusion_baseline"
)

CHECKPOINT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

RESULT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


def set_seed(seed=SEED):

    random.seed(seed)
    np.random.seed(seed)

    torch.manual_seed(seed)

    if torch.cuda.is_available():
        torch.cuda.manual_seed_all(seed)


def load_features(split):

    path = FEATURE_ROOT / f"{split}.pt"

    data = torch.load(
        path,
        map_location="cpu",
        weights_only=False
    )

    return data


def standardize(
    train,
    validation,
    test
):

    mean = train.mean(
        dim=0,
        keepdim=True
    )

    std = train.std(
        dim=0,
        keepdim=True
    )

    std = torch.where(
        std < 1e-6,
        torch.ones_like(std),
        std
    )

    train = (
        train - mean
    ) / std

    validation = (
        validation - mean
    ) / std

    test = (
        test - mean
    ) / std

    return (
        train,
        validation,
        test,
        mean,
        std
    )


class FusionMLP(nn.Module):

    def __init__(
        self,
        input_dim=2816
    ):

        super().__init__()

        self.network = nn.Sequential(

            nn.Linear(
                input_dim,
                512
            ),

            nn.ReLU(),

            nn.Dropout(
                0.30
            ),

            nn.Linear(
                512,
                128
            ),

            nn.ReLU(),

            nn.Dropout(
                0.20
            ),

            nn.Linear(
                128,
                2
            )
        )

    def forward(self, x):

        return self.network(x)


# END REGISTERED SOURCE BLOCK


In [26]:
%%project_source multimodal-fake-news-detection/scripts/train_multimodal_fusion.py 1
def compute_metrics(
    labels,
    predictions,
    probabilities
):

    metrics = {

        "accuracy":
            accuracy_score(
                labels,
                predictions
            ),

        "precision":
            precision_score(
                labels,
                predictions,
                zero_division=0
            ),

        "recall":
            recall_score(
                labels,
                predictions,
                zero_division=0
            ),

        "f1":
            f1_score(
                labels,
                predictions,
                zero_division=0
            ),

        "f1_macro":
            f1_score(
                labels,
                predictions,
                average="macro",
                zero_division=0
            ),
    }

    try:

        metrics["roc_auc"] = (
            roc_auc_score(
                labels,
                probabilities
            )
        )

    except ValueError:

        metrics["roc_auc"] = None


    try:

        metrics["pr_auc"] = (
            average_precision_score(
                labels,
                probabilities
            )
        )

    except ValueError:

        metrics["pr_auc"] = None


    return metrics


def evaluate(
    model,
    loader,
    criterion,
    device
):

    model.eval()

    total_loss = 0.0

    labels_all = []
    predictions_all = []
    probabilities_all = []

    with torch.no_grad():

        for features, labels in loader:

            features = features.to(
                device,
                non_blocking=True
            )

            labels = labels.to(
                device,
                non_blocking=True
            )

            logits = model(
                features
            )

            loss = criterion(
                logits,
                labels
            )

            probabilities = (
                torch.softmax(
                    logits,
                    dim=1
                )[:, 1]
            )

            predictions = (
                torch.argmax(
                    logits,
                    dim=1
                )
            )

            total_loss += (
                loss.item()
            )

            labels_all.extend(
                labels.cpu()
                .numpy()
                .tolist()
            )

            predictions_all.extend(
                predictions.cpu()
                .numpy()
                .tolist()
            )

            probabilities_all.extend(
                probabilities.cpu()
                .numpy()
                .tolist()
            )


    metrics = compute_metrics(
        labels_all,
        predictions_all,
        probabilities_all
    )

    metrics["loss"] = (
        total_loss
        / len(loader)
    )

    return (
        metrics,
        labels_all,
        predictions_all,
        probabilities_all
    )


# END REGISTERED SOURCE BLOCK


In [27]:
%%project_source multimodal-fake-news-detection/scripts/train_multimodal_fusion.py 2
def train_epoch(
    model,
    loader,
    optimizer,
    criterion,
    device
):

    model.train()

    total_loss = 0.0

    for features, labels in loader:

        features = features.to(
            device,
            non_blocking=True
        )

        labels = labels.to(
            device,
            non_blocking=True
        )

        optimizer.zero_grad(
            set_to_none=True
        )

        logits = model(
            features
        )

        loss = criterion(
            logits,
            labels
        )

        loss.backward()

        torch.nn.utils.clip_grad_norm_(
            model.parameters(),
            max_norm=1.0
        )

        optimizer.step()

        total_loss += (
            loss.item()
        )

    return (
        total_loss / len(loader)
    )


def main():

    parser = argparse.ArgumentParser()

    parser.add_argument(
        "--epochs",
        type=int,
        default=30
    )

    parser.add_argument(
        "--batch-size",
        type=int,
        default=256
    )

    parser.add_argument(
        "--lr",
        type=float,
        default=1e-3
    )

    parser.add_argument(
        "--smoke-test",
        action="store_true"
    )

    args = parser.parse_args()

    set_seed()

    device = torch.device(
        "cuda"
        if torch.cuda.is_available()
        else "cpu"
    )


    print("=" * 70)
    print("MULTIMODAL FUSION BASELINE")
    print("=" * 70)

    print(
        f"\nDevice: {device}"
    )

    if device.type == "cuda":

        print(
            "GPU:",
            torch.cuda.get_device_name(0)
        )


    # --------------------------------------------------------
    # Load extracted features
    # --------------------------------------------------------

    train = load_features(
        "train"
    )

    validation = load_features(
        "validation"
    )

    test = load_features(
        "test"
    )


    train_text = (
        train["text_features"]
        .float()
    )

    validation_text = (
        validation["text_features"]
        .float()
    )

    test_text = (
        test["text_features"]
        .float()
    )


    train_image = (
        train["image_features"]
        .float()
    )

    validation_image = (
        validation["image_features"]
        .float()
    )

    test_image = (
        test["image_features"]
        .float()
    )


    # --------------------------------------------------------
    # Normalize each modality independently.
    # Statistics are estimated from TRAIN ONLY.
    # --------------------------------------------------------

    (
        train_text,
        validation_text,
        test_text,
        text_mean,
        text_std
    ) = standardize(
        train_text,
        validation_text,
        test_text
    )


    (
        train_image,
        validation_image,
        test_image,
        image_mean,
        image_std
    ) = standardize(
        train_image,
        validation_image,
        test_image
    )


    # --------------------------------------------------------
    # Concatenate modalities
    # --------------------------------------------------------

    train_features = torch.cat(
        [
            train_text,
            train_image
        ],
        dim=1
    )

    validation_features = torch.cat(
        [
            validation_text,
            validation_image
        ],
        dim=1
    )

    test_features = torch.cat(
        [
            test_text,
            test_image
        ],
        dim=1
    )


    train_labels = (
        train["labels"].long()
    )

    validation_labels = (
        validation["labels"].long()
    )

    test_labels = (
        test["labels"].long()
    )


    train_ids = train["ids"]
    validation_ids = validation["ids"]
    test_ids = test["ids"]


    print("\nFeature shapes:")

    print(
        "Train:     ",
        tuple(
            train_features.shape
        )
    )

    print(
        "Validation:",
        tuple(
            validation_features.shape
        )
    )

    print(
        "Test:      ",
        tuple(
            test_features.shape
        )
    )


    if (
        train_features.shape[1]
        != 2816
    ):

        raise ValueError(
            "Expected 2816 fused features."
        )


    # --------------------------------------------------------
    # Smoke test
    # --------------------------------------------------------

    if args.smoke_test:

        print(
            "\nSMOKE TEST MODE"
        )

        train_features = (
            train_features[:512]
        )

        train_labels = (
            train_labels[:512]
        )

        train_ids = (
            train_ids[:512]
        )

        validation_features = (
            validation_features[:256]
        )

        validation_labels = (
            validation_labels[:256]
        )

        validation_ids = (
            validation_ids[:256]
        )

        test_features = (
            test_features[:256]
        )

        test_labels = (
            test_labels[:256]
        )

        test_ids = (
            test_ids[:256]
        )

        args.epochs = 3


    print("\nDataset sizes:")

    print(
        f"Train:      "
        f"{len(train_labels):,}"
    )

    print(
        f"Validation: "
        f"{len(validation_labels):,}"
    )

    print(
        f"Test:       "
        f"{len(test_labels):,}"
    )


    train_dataset = TensorDataset(
        train_features,
        train_labels
    )

    validation_dataset = TensorDataset(
        validation_features,
        validation_labels
    )

    test_dataset = TensorDataset(
        test_features,
        test_labels
    )


    train_loader = DataLoader(
        train_dataset,
        batch_size=args.batch_size,
        shuffle=True,
        pin_memory=(
            device.type == "cuda"
        )
    )

    validation_loader = DataLoader(
        validation_dataset,
        batch_size=args.batch_size,
        shuffle=False,
        pin_memory=(
            device.type == "cuda"
        )
    )

    test_loader = DataLoader(
        test_dataset,
        batch_size=args.batch_size,
        shuffle=False,
        pin_memory=(
            device.type == "cuda"
        )
    )


    model = FusionMLP().to(
        device
    )


    criterion = (
        nn.CrossEntropyLoss()
    )


    optimizer = AdamW(
        model.parameters(),
        lr=args.lr,
        weight_decay=1e-4
    )


    best_macro_f1 = -1.0
    epochs_without_improvement = 0
    patience = 5

    history = []


    # --------------------------------------------------------
    # Training
    # --------------------------------------------------------

    for epoch in range(
        1,
        args.epochs + 1
    ):

        print(
            "\n" + "=" * 70
        )

        print(
            f"EPOCH "
            f"{epoch}/{args.epochs}"
        )

        print("=" * 70)


        train_loss = train_epoch(
            model,
            train_loader,
            optimizer,
            criterion,
            device
        )


        (
            validation_metrics,
            _,
            _,
            _
        ) = evaluate(
            model,
            validation_loader,
            criterion,
            device
        )


        print(
            f"\nTrain loss: "
            f"{train_loss:.4f}"
        )


        print(
            "\nValidation metrics:"
        )


        for name, value in (
            validation_metrics.items()
        ):

            if value is None:

                print(
                    f"{name:12s}: N/A"
                )

            else:

                print(
                    f"{name:12s}: "
                    f"{value:.4f}"
                )


        history.append({

            "epoch":
                epoch,

            "train_loss":
                train_loss,

            **{
                f"validation_{k}":
                    v

                for k, v
                in validation_metrics.items()
            }
        })


        current_macro_f1 = (
            validation_metrics[
                "f1_macro"
            ]
        )


        if (
            current_macro_f1
            > best_macro_f1
        ):

            best_macro_f1 = (
                current_macro_f1
            )

            epochs_without_improvement = 0

            print(
                "\nNew best validation "
                "macro F1. "
                "Saving checkpoint."
            )


            torch.save(
                {
                    "model_state_dict":
                        model.state_dict(),

                    "text_mean":
                        text_mean,

                    "text_std":
                        text_std,

                    "image_mean":
                        image_mean,

                    "image_std":
                        image_std,

                    "validation_macro_f1":
                        best_macro_f1,

                    "input_dim":
                        2816,
                },

                CHECKPOINT_ROOT
                / "best_model.pt"
            )


        else:

            epochs_without_improvement += 1

            print(
                "\nNo validation macro "
                "F1 improvement."
            )


            if (
                epochs_without_improvement
                >= patience
            ):

                print(
                    "Early stopping "
                    "triggered."
                )

                break


    # --------------------------------------------------------
    # Save history
    # --------------------------------------------------------

    pd.DataFrame(
        history
    ).to_csv(
        RESULT_ROOT
        / "training_history.csv",
        index=False
    )


    # --------------------------------------------------------
    # Load best fusion model
    # --------------------------------------------------------

    print(
        "\nLoading best checkpoint..."
    )


    checkpoint = torch.load(
        CHECKPOINT_ROOT
        / "best_model.pt",
        map_location=device,
        weights_only=False
    )


    model.load_state_dict(
        checkpoint[
            "model_state_dict"
        ]
    )


    # --------------------------------------------------------
    # Test evaluation
    # --------------------------------------------------------

    (
        test_metrics,
        labels,
        predictions,
        probabilities
    ) = evaluate(
        model,
        test_loader,
        criterion,
        device
    )


    print(
        "\n" + "=" * 70
    )

    print(
        "TEST RESULTS"
    )

    print("=" * 70)


    for name, value in (
        test_metrics.items()
    ):

        if value is None:

            print(
                f"{name:12s}: N/A"
            )

        else:

            print(
                f"{name:12s}: "
                f"{value:.4f}"
            )


    matrix = confusion_matrix(
        labels,
        predictions
    )


    print(
        "\nConfusion matrix:"
    )

    print(matrix)


    # --------------------------------------------------------
    # Save results
    # --------------------------------------------------------

    with (
        RESULT_ROOT
        / "test_metrics.json"
    ).open(
        "w",
        encoding="utf-8"
    ) as f:

        json.dump(
            {
                **test_metrics,

                "confusion_matrix":
                    matrix.tolist(),

                "best_validation_macro_f1":
                    best_macro_f1,

                "model":
                    "frozen_feature_concat_mlp",

                "text_encoder":
                    "fine_tuned_roberta_base",

                "image_encoder":
                    "fine_tuned_resnet50",

                "text_dimension":
                    768,

                "image_dimension":
                    2048,

                "fusion_dimension":
                    2816,

                "seed":
                    SEED,

                "batch_size":
                    args.batch_size,

                "learning_rate":
                    args.lr,
            },

            f,
            indent=2
        )


    prediction_df = pd.DataFrame({

        "id":
            test_ids,

        "label":
            labels,

        "prediction":
            predictions,

        "probability_class_1":
            probabilities
    })


    prediction_df.to_csv(
        RESULT_ROOT
        / "test_predictions.csv",
        index=False
    )


    print(
        "\nResults saved to:",
        RESULT_ROOT
    )

    print(
        "Best model saved to:",
        CHECKPOINT_ROOT
    )


# END REGISTERED SOURCE BLOCK


In [28]:
%%project_source multimodal-fake-news-detection/scripts/train_multimodal_fusion.py 3
if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


### 5.3 Tune multimodal fusion

Compare development fusion settings to investigate generalisation and overfitting; these are development experiments.

**Source:** `multimodal-fake-news-detection/scripts/tune_multimodal_fusion.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `random`, `sklearn`, `torch`  
**Top-level components:** `set_seed`, `load_split`, `standardise`, `FusionMLP`, `evaluate`, `run_experiment`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/multimodal_features`
- `results/metrics/multimodal_fusion_tuning`

The following cells contain the complete source; Run All registers it for inspection/export.

In [29]:
%%project_source multimodal-fake-news-detection/scripts/tune_multimodal_fusion.py 0
import json
import random
from pathlib import Path

import numpy as np
import pandas as pd
import torch
import torch.nn as nn

from torch.utils.data import (
    DataLoader,
    TensorDataset,
)

from sklearn.metrics import (
    accuracy_score,
    f1_score,
)


FEATURE_ROOT = Path(
    "data/processed/fakeddit/multimodal_features"
)

OUTPUT_ROOT = Path(
    "results/metrics/multimodal_fusion_tuning"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


SEEDS = [42, 52, 62]

MAX_EPOCHS = 25
PATIENCE = 4
BATCH_SIZE = 256


CONFIGS = [
    {
        "name": "bottleneck_64",
        "hidden": [64],
        "dropout": [0.30],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        "name": "small_128",
        "hidden": [128],
        "dropout": [0.30],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        "name": "small_128_high_dropout",
        "hidden": [128],
        "dropout": [0.50],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        "name": "medium_256",
        "hidden": [256],
        "dropout": [0.30],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        "name": "medium_256_high_dropout",
        "hidden": [256],
        "dropout": [0.50],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        "name": "two_layer_128_64",
        "hidden": [128, 64],
        "dropout": [0.40, 0.30],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        "name": "two_layer_256_64",
        "hidden": [256, 64],
        "dropout": [0.40, 0.30],
        "lr": 3e-4,
        "weight_decay": 1e-3,
    },

    {
        # Similar to the previous high-capacity baseline,
        # included as a control.
        "name": "large_512_128",
        "hidden": [512, 128],
        "dropout": [0.30, 0.20],
        "lr": 1e-3,
        "weight_decay": 1e-4,
    },
]


def set_seed(seed):

    random.seed(seed)
    np.random.seed(seed)

    torch.manual_seed(seed)

    if torch.cuda.is_available():

        torch.cuda.manual_seed_all(
            seed
        )


def load_split(split):

    data = torch.load(
        FEATURE_ROOT / f"{split}.pt",
        map_location="cpu",
        weights_only=False
    )

    text = (
        data["text_features"]
        .float()
    )

    image = (
        data["image_features"]
        .float()
    )

    labels = (
        data["labels"]
        .long()
    )

    return (
        text,
        image,
        labels
    )


def standardise(
    train_tensor,
    validation_tensor
):

    mean = train_tensor.mean(
        dim=0,
        keepdim=True
    )

    std = train_tensor.std(
        dim=0,
        keepdim=True
    )

    std = torch.where(
        std < 1e-6,
        torch.ones_like(std),
        std
    )

    train_scaled = (
        train_tensor - mean
    ) / std

    validation_scaled = (
        validation_tensor - mean
    ) / std

    return (
        train_scaled,
        validation_scaled
    )


# END REGISTERED SOURCE BLOCK


In [30]:
%%project_source multimodal-fake-news-detection/scripts/tune_multimodal_fusion.py 1
class FusionMLP(nn.Module):

    def __init__(
        self,
        input_dim,
        hidden_dims,
        dropout_values
    ):

        super().__init__()

        layers = []

        current_dim = input_dim

        for hidden_dim, dropout in zip(
            hidden_dims,
            dropout_values
        ):

            layers.extend([
                nn.Linear(
                    current_dim,
                    hidden_dim
                ),

                nn.ReLU(),

                nn.Dropout(
                    dropout
                ),
            ])

            current_dim = hidden_dim

        layers.append(
            nn.Linear(
                current_dim,
                2
            )
        )

        self.network = nn.Sequential(
            *layers
        )

    def forward(self, x):

        return self.network(x)


@torch.no_grad()
def evaluate(
    model,
    loader,
    criterion,
    device
):

    model.eval()

    losses = []

    labels_all = []
    predictions_all = []

    for features, labels in loader:

        features = features.to(
            device,
            non_blocking=True
        )

        labels = labels.to(
            device,
            non_blocking=True
        )

        logits = model(
            features
        )

        loss = criterion(
            logits,
            labels
        )

        losses.append(
            loss.item()
            * labels.size(0)
        )

        predictions = torch.argmax(
            logits,
            dim=1
        )

        labels_all.extend(
            labels.cpu().numpy()
        )

        predictions_all.extend(
            predictions.cpu().numpy()
        )

    labels_all = np.asarray(
        labels_all
    )

    predictions_all = np.asarray(
        predictions_all
    )

    return {
        "loss":
            float(
                sum(losses)
                / len(labels_all)
            ),

        "accuracy":
            float(
                accuracy_score(
                    labels_all,
                    predictions_all
                )
            ),

        "f1_macro":
            float(
                f1_score(
                    labels_all,
                    predictions_all,
                    average="macro"
                )
            ),
    }


def run_experiment(
    config,
    seed,
    train_loader,
    validation_loader,
    input_dim,
    device
):

    set_seed(seed)

    model = FusionMLP(
        input_dim=input_dim,
        hidden_dims=config["hidden"],
        dropout_values=config["dropout"]
    ).to(device)

    criterion = (
        nn.CrossEntropyLoss()
    )

    optimizer = torch.optim.AdamW(
        model.parameters(),
        lr=config["lr"],
        weight_decay=config[
            "weight_decay"
        ]
    )

    best_macro_f1 = -1.0
    best_epoch = None
    best_accuracy = None
    best_loss = None

    epochs_without_improvement = 0

    for epoch in range(
        1,
        MAX_EPOCHS + 1
    ):

        model.train()

        for features, labels in train_loader:

            features = features.to(
                device,
                non_blocking=True
            )

            labels = labels.to(
                device,
                non_blocking=True
            )

            optimizer.zero_grad(
                set_to_none=True
            )

            logits = model(
                features
            )

            loss = criterion(
                logits,
                labels
            )

            loss.backward()

            torch.nn.utils.clip_grad_norm_(
                model.parameters(),
                max_norm=1.0
            )

            optimizer.step()

        validation_metrics = evaluate(
            model,
            validation_loader,
            criterion,
            device
        )

        macro_f1 = (
            validation_metrics[
                "f1_macro"
            ]
        )

        if (
            macro_f1
            > best_macro_f1 + 1e-5
        ):

            best_macro_f1 = (
                macro_f1
            )

            best_epoch = epoch

            best_accuracy = (
                validation_metrics[
                    "accuracy"
                ]
            )

            best_loss = (
                validation_metrics[
                    "loss"
                ]
            )

            epochs_without_improvement = 0

        else:

            epochs_without_improvement += 1

        if (
            epochs_without_improvement
            >= PATIENCE
        ):
            break

    return {
        "config":
            config["name"],

        "seed":
            seed,

        "best_epoch":
            int(best_epoch),

        "validation_macro_f1":
            float(best_macro_f1),

        "validation_accuracy":
            float(best_accuracy),

        "validation_loss":
            float(best_loss),
    }


# END REGISTERED SOURCE BLOCK


In [31]:
%%project_source multimodal-fake-news-detection/scripts/tune_multimodal_fusion.py 2
def main():

    device = torch.device(
        "cuda"
        if torch.cuda.is_available()
        else "cpu"
    )

    print("=" * 70)
    print("MULTIMODAL FUSION TUNING")
    print("=" * 70)

    print(
        f"\nDevice: {device}"
    )

    if device.type == "cuda":

        print(
            "GPU:",
            torch.cuda.get_device_name(0)
        )


    # --------------------------------------------------------
    # TRAIN + VALIDATION ONLY
    # --------------------------------------------------------

    train_text, train_image, train_labels = (
        load_split("train")
    )

    validation_text, validation_image, validation_labels = (
        load_split("validation")
    )


    # Standardise each modality separately.
    # Statistics are learned from TRAIN only.
    train_text, validation_text = (
        standardise(
            train_text,
            validation_text
        )
    )

    train_image, validation_image = (
        standardise(
            train_image,
            validation_image
        )
    )


    train_features = torch.cat(
        [
            train_text,
            train_image
        ],
        dim=1
    )

    validation_features = torch.cat(
        [
            validation_text,
            validation_image
        ],
        dim=1
    )


    print(
        "\nTraining samples:",
        len(train_labels)
    )

    print(
        "Validation samples:",
        len(validation_labels)
    )

    print(
        "Feature dimension:",
        train_features.shape[1]
    )

    print(
        "\nTEST SET IS NOT LOADED."
    )


    train_dataset = TensorDataset(
        train_features,
        train_labels
    )

    validation_dataset = TensorDataset(
        validation_features,
        validation_labels
    )


    validation_loader = DataLoader(
        validation_dataset,
        batch_size=BATCH_SIZE,
        shuffle=False,
        pin_memory=(
            device.type == "cuda"
        )
    )


    all_runs = []


    for config in CONFIGS:

        print(
            "\n" + "=" * 70
        )

        print(
            config["name"].upper()
        )

        print("=" * 70)

        print(
            "Hidden:",
            config["hidden"]
        )

        print(
            "Dropout:",
            config["dropout"]
        )

        print(
            "LR:",
            config["lr"]
        )

        print(
            "Weight decay:",
            config["weight_decay"]
        )


        for seed in SEEDS:

            # Recreate shuffled loader
            # using this experiment's seed.
            generator = (
                torch.Generator()
            )

            generator.manual_seed(
                seed
            )

            train_loader = DataLoader(
                train_dataset,
                batch_size=BATCH_SIZE,
                shuffle=True,
                generator=generator,
                pin_memory=(
                    device.type == "cuda"
                )
            )


            result = run_experiment(
                config=config,
                seed=seed,
                train_loader=train_loader,
                validation_loader=validation_loader,
                input_dim=(
                    train_features.shape[1]
                ),
                device=device
            )

            all_runs.append(
                result
            )

            print(
                f"Seed {seed}: "
                f"best epoch "
                f"{result['best_epoch']:2d} | "
                f"macro F1 "
                f"{result['validation_macro_f1']:.4f} | "
                f"accuracy "
                f"{result['validation_accuracy']:.4f}"
            )


    runs_df = pd.DataFrame(
        all_runs
    )

    runs_df.to_csv(
        OUTPUT_ROOT
        / "all_runs.csv",
        index=False
    )


    summary = (
        runs_df
        .groupby("config")
        .agg(
            mean_macro_f1=(
                "validation_macro_f1",
                "mean"
            ),

            std_macro_f1=(
                "validation_macro_f1",
                "std"
            ),

            mean_accuracy=(
                "validation_accuracy",
                "mean"
            ),

            mean_best_epoch=(
                "best_epoch",
                "mean"
            ),
        )
        .sort_values(
            "mean_macro_f1",
            ascending=False
        )
        .reset_index()
    )


    summary.to_csv(
        OUTPUT_ROOT
        / "summary.csv",
        index=False
    )


    print(
        "\n" + "=" * 70
    )

    print(
        "VALIDATION-ONLY RANKING"
    )

    print("=" * 70)

    print(
        summary.to_string(
            index=False,
            float_format=lambda x:
                f"{x:.4f}"
        )
    )


    best_name = (
        summary.iloc[0][
            "config"
        ]
    )

    best_config = next(
        config
        for config in CONFIGS
        if config["name"]
        == best_name
    )


    best_result = {
        "selection_metric":
            "mean validation macro F1",

        "seeds":
            SEEDS,

        "test_evaluated":
            False,

        "best_config":
            best_config,

        "validation_summary":
            summary.iloc[0]
            .to_dict(),
    }


    with (
        OUTPUT_ROOT
        / "best_config.json"
    ).open(
        "w",
        encoding="utf-8"
    ) as f:

        json.dump(
            best_result,
            f,
            indent=2
        )


    print(
        "\nSelected configuration:"
    )

    print(
        json.dumps(
            best_config,
            indent=2
        )
    )

    print(
        "\nNo test evaluation "
        "was performed."
    )

    print(
        "\nResults saved to:",
        OUTPUT_ROOT
    )


# END REGISTERED SOURCE BLOCK


In [32]:
%%project_source multimodal-fake-news-detection/scripts/tune_multimodal_fusion.py 3
if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


### 5.4 Evaluate linear fusion

Compare linear probes over text, image and combined representations as a simpler fusion control.

**Source:** `multimodal-fake-news-detection/scripts/evaluate_linear_fusion.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `sklearn`, `torch`  
**Top-level components:** `load_split`, `metrics`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/multimodal_features`
- `results/metrics/linear_fusion_ablation`

The following cells contain the complete source; Run All registers it for inspection/export.

In [33]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_linear_fusion.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd
import torch

from sklearn.linear_model import LogisticRegression
from sklearn.preprocessing import StandardScaler
from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
    confusion_matrix,
)


FEATURE_ROOT = Path(
    "data/processed/fakeddit/multimodal_features"
)

RESULT_ROOT = Path(
    "results/metrics/linear_fusion_ablation"
)

RESULT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

SEED = 42


def load_split(split):

    data = torch.load(
        FEATURE_ROOT / f"{split}.pt",
        map_location="cpu",
        weights_only=False
    )

    return {
        "ids": list(data["ids"]),
        "labels": data["labels"].numpy(),
        "text": data["text_features"].numpy(),
        "image": data["image_features"].numpy(),
    }


def metrics(
    y_true,
    y_pred,
    y_prob
):

    return {
        "accuracy": float(
            accuracy_score(
                y_true,
                y_pred
            )
        ),

        "precision": float(
            precision_score(
                y_true,
                y_pred,
                zero_division=0
            )
        ),

        "recall": float(
            recall_score(
                y_true,
                y_pred,
                zero_division=0
            )
        ),

        "f1": float(
            f1_score(
                y_true,
                y_pred,
                zero_division=0
            )
        ),

        "f1_macro": float(
            f1_score(
                y_true,
                y_pred,
                average="macro",
                zero_division=0
            )
        ),

        "roc_auc": float(
            roc_auc_score(
                y_true,
                y_prob
            )
        ),

        "pr_auc": float(
            average_precision_score(
                y_true,
                y_prob
            )
        ),

        "confusion_matrix":
            confusion_matrix(
                y_true,
                y_pred
            ).tolist(),
    }


train = load_split("train")
validation = load_split("validation")
test = load_split("test")


experiments = {
    "text_only": (
        train["text"],
        validation["text"],
        test["text"]
    ),

    "image_only": (
        train["image"],
        validation["image"],
        test["image"]
    ),

    "text_image_concat": (
        np.concatenate(
            [
                train["text"],
                train["image"]
            ],
            axis=1
        ),

        np.concatenate(
            [
                validation["text"],
                validation["image"]
            ],
            axis=1
        ),

        np.concatenate(
            [
                test["text"],
                test["image"]
            ],
            axis=1
        ),
    )
}


# END REGISTERED SOURCE BLOCK


In [34]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_linear_fusion.py 1
all_results = {}


for name, (
    X_train,
    X_validation,
    X_test
) in experiments.items():

    print("\n" + "=" * 70)
    print(name.upper())
    print("=" * 70)

    print(
        "Dimensions:",
        X_train.shape[1]
    )

    # Fit scaling using TRAIN ONLY.
    scaler = StandardScaler()

    X_train = scaler.fit_transform(
        X_train
    )

    X_validation = scaler.transform(
        X_validation
    )

    X_test = scaler.transform(
        X_test
    )


    model = LogisticRegression(
        C=1.0,
        max_iter=3000,
        solver="lbfgs",
        random_state=SEED
    )


    print("Training...")

    model.fit(
        X_train,
        train["labels"]
    )


    # --------------------------------------------------------
    # Validation
    # --------------------------------------------------------

    validation_prob = (
        model.predict_proba(
            X_validation
        )[:, 1]
    )

    validation_pred = (
        model.predict(
            X_validation
        )
    )

    validation_metrics = metrics(
        validation["labels"],
        validation_pred,
        validation_prob
    )


    print(
        "\nValidation metrics:"
    )

    for key, value in (
        validation_metrics.items()
    ):

        if key == "confusion_matrix":
            continue

        print(
            f"{key:12s}: "
            f"{value:.4f}"
        )


    print(
        "Confusion matrix:"
    )

    print(
        np.array(
            validation_metrics[
                "confusion_matrix"
            ]
        )
    )


    # --------------------------------------------------------
    # Test
    # --------------------------------------------------------

    test_prob = (
        model.predict_proba(
            X_test
        )[:, 1]
    )

    test_pred = (
        model.predict(
            X_test
        )
    )

    test_metrics = metrics(
        test["labels"],
        test_pred,
        test_prob
    )


    print(
        "\nTest metrics:"
    )

    for key, value in (
        test_metrics.items()
    ):

        if key == "confusion_matrix":
            continue

        print(
            f"{key:12s}: "
            f"{value:.4f}"
        )


    print(
        "Confusion matrix:"
    )

    print(
        np.array(
            test_metrics[
                "confusion_matrix"
            ]
        )
    )


    all_results[name] = {
        "validation":
            validation_metrics,

        "test":
            test_metrics,

        "feature_dimension":
            int(X_train.shape[1]),

        "classifier":
            "logistic_regression",

        "C":
            1.0
    }


    predictions = pd.DataFrame({
        "id":
            test["ids"],

        "label":
            test["labels"],

        "prediction":
            test_pred,

        "probability_class_1":
            test_prob
    })


    predictions.to_csv(
        RESULT_ROOT
        / f"{name}_test_predictions.csv",
        index=False
    )


# END REGISTERED SOURCE BLOCK


In [35]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_linear_fusion.py 2
with (
    RESULT_ROOT
    / "results.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        all_results,
        f,
        indent=2
    )


print("\n" + "=" * 70)
print("LINEAR FUSION ABLATION COMPLETE")
print("=" * 70)

print(
    "\nResults saved to:",
    RESULT_ROOT
)
# END REGISTERED SOURCE BLOCK


### 5.5 Export baseline probabilities

Run the locked unimodal checkpoints and export per-ID class probabilities for paired fusion.

**Source:** `multimodal-fake-news-detection/scripts/export_baseline_probabilities.py`  
**Imported modules:** `PIL`, `pandas`, `pathlib`, `torch`, `torchvision`, `transformers`  
**Top-level components:** `TextDataset`, `ImageDataset`, `export_roberta`, `export_resnet`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/development_clean`
- `checkpoints/roberta_baseline`
- `checkpoints/resnet50_baseline/best_model.pt`
- `results/metrics/baseline_probabilities`

The following cells contain the complete source; Run All registers it for inspection/export.

In [36]:
%%project_source multimodal-fake-news-detection/scripts/export_baseline_probabilities.py 0
from pathlib import Path

import pandas as pd
from PIL import Image

import torch
import torch.nn as nn
from torch.utils.data import Dataset, DataLoader

from transformers import (
    AutoTokenizer,
    AutoModelForSequenceClassification,
)

from torchvision.models import resnet50
from torchvision import transforms


DATA_ROOT = Path(
    "data/processed/fakeddit/development_clean"
)

ROBERTA_CHECKPOINT = Path(
    "checkpoints/roberta_baseline"
)

RESNET_CHECKPOINT = Path(
    "checkpoints/resnet50_baseline/best_model.pt"
)

OUTPUT_ROOT = Path(
    "results/metrics/baseline_probabilities"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

MAX_LENGTH = 64
BATCH_SIZE_TEXT = 16
BATCH_SIZE_IMAGE = 32
NUM_WORKERS = 4


class TextDataset(Dataset):

    def __init__(
        self,
        dataframe,
        tokenizer
    ):

        self.df = (
            dataframe
            .reset_index(drop=True)
        )

        self.tokenizer = tokenizer

    def __len__(self):
        return len(self.df)

    def __getitem__(self, idx):

        row = self.df.iloc[idx]

        tokens = self.tokenizer(
            str(row["text"]),
            padding="max_length",
            truncation=True,
            max_length=MAX_LENGTH,
            return_tensors="pt"
        )

        return {
            "id": str(row["id"]),

            "label": int(
                row["label"]
            ),

            "input_ids":
                tokens["input_ids"]
                .squeeze(0),

            "attention_mask":
                tokens["attention_mask"]
                .squeeze(0),
        }


class ImageDataset(Dataset):

    def __init__(
        self,
        dataframe,
        transform
    ):

        self.df = (
            dataframe
            .reset_index(drop=True)
        )

        self.transform = transform

    def __len__(self):
        return len(self.df)

    def __getitem__(self, idx):

        row = self.df.iloc[idx]

        image_path = Path(
            str(row["image_path"])
        )

        with Image.open(
            image_path
        ) as image:

            image = image.convert(
                "RGB"
            )

            image = self.transform(
                image
            )

        return {
            "id": str(row["id"]),

            "label": int(
                row["label"]
            ),

            "image": image,
        }


@torch.no_grad()
def export_roberta(
    dataframe,
    split,
    model,
    tokenizer,
    device
):

    dataset = TextDataset(
        dataframe,
        tokenizer
    )

    loader = DataLoader(
        dataset,
        batch_size=BATCH_SIZE_TEXT,
        shuffle=False,
        num_workers=0,
        pin_memory=(
            device.type == "cuda"
        )
    )

    ids = []
    labels = []
    probabilities = []
    predictions = []

    model.eval()

    for batch in loader:

        input_ids = (
            batch["input_ids"]
            .to(
                device,
                non_blocking=True
            )
        )

        attention_mask = (
            batch["attention_mask"]
            .to(
                device,
                non_blocking=True
            )
        )

        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=(
                device.type == "cuda"
            )
        ):

            outputs = model(
                input_ids=input_ids,
                attention_mask=attention_mask
            )

            logits = outputs.logits

        probs = torch.softmax(
            logits,
            dim=1
        )[:, 1]

        preds = torch.argmax(
            logits,
            dim=1
        )

        ids.extend(
            batch["id"]
        )

        labels.extend(
            batch["label"]
            .numpy()
            .tolist()
        )

        probabilities.extend(
            probs
            .cpu()
            .numpy()
            .tolist()
        )

        predictions.extend(
            preds
            .cpu()
            .numpy()
            .tolist()
        )

    output = pd.DataFrame({
        "id": ids,
        "label": labels,
        "prediction": predictions,
        "probability_class_1":
            probabilities,
    })

    path = (
        OUTPUT_ROOT
        / f"roberta_{split}.csv"
    )

    output.to_csv(
        path,
        index=False
    )

    print(
        f"RoBERTa {split}: "
        f"{len(output):,} rows -> {path}"
    )


# END REGISTERED SOURCE BLOCK


In [37]:
%%project_source multimodal-fake-news-detection/scripts/export_baseline_probabilities.py 1
@torch.no_grad()
def export_resnet(
    dataframe,
    split,
    model,
    transform,
    device
):

    dataset = ImageDataset(
        dataframe,
        transform
    )

    loader_kwargs = {
        "batch_size":
            BATCH_SIZE_IMAGE,

        "shuffle":
            False,

        "num_workers":
            NUM_WORKERS,

        "pin_memory":
            device.type == "cuda",
    }

    if NUM_WORKERS > 0:
        loader_kwargs[
            "persistent_workers"
        ] = True

    loader = DataLoader(
        dataset,
        **loader_kwargs
    )

    ids = []
    labels = []
    probabilities = []
    predictions = []

    model.eval()

    for batch in loader:

        images = (
            batch["image"]
            .to(
                device,
                non_blocking=True
            )
        )

        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=(
                device.type == "cuda"
            )
        ):

            logits = model(
                images
            )

        probs = torch.softmax(
            logits,
            dim=1
        )[:, 1]

        preds = torch.argmax(
            logits,
            dim=1
        )

        ids.extend(
            batch["id"]
        )

        labels.extend(
            batch["label"]
            .numpy()
            .tolist()
        )

        probabilities.extend(
            probs
            .cpu()
            .numpy()
            .tolist()
        )

        predictions.extend(
            preds
            .cpu()
            .numpy()
            .tolist()
        )

    output = pd.DataFrame({
        "id": ids,
        "label": labels,
        "prediction": predictions,
        "probability_class_1":
            probabilities,
    })

    path = (
        OUTPUT_ROOT
        / f"resnet_{split}.csv"
    )

    output.to_csv(
        path,
        index=False
    )

    print(
        f"ResNet {split}: "
        f"{len(output):,} rows -> {path}"
    )


def main():

    device = torch.device(
        "cuda"
        if torch.cuda.is_available()
        else "cpu"
    )

    print("=" * 70)
    print("EXPORT BASELINE PROBABILITIES")
    print("=" * 70)

    print(
        f"\nDevice: {device}"
    )

    if device.type == "cuda":

        print(
            "GPU:",
            torch.cuda.get_device_name(0)
        )


    # --------------------------------------------------------
    # RoBERTa
    # --------------------------------------------------------

    print(
        "\nLoading RoBERTa checkpoint..."
    )

    tokenizer = (
        AutoTokenizer
        .from_pretrained(
            ROBERTA_CHECKPOINT
        )
    )

    roberta = (
        AutoModelForSequenceClassification
        .from_pretrained(
            ROBERTA_CHECKPOINT
        )
    )

    roberta.to(device)


    # --------------------------------------------------------
    # ResNet
    # --------------------------------------------------------

    print(
        "Loading ResNet checkpoint..."
    )

    resnet_checkpoint = torch.load(
        RESNET_CHECKPOINT,
        map_location="cpu",
        weights_only=True
    )

    resnet = resnet50(
        weights=None
    )

    features = (
        resnet.fc.in_features
    )

    resnet.fc = nn.Linear(
        features,
        2
    )

    resnet.load_state_dict(
        resnet_checkpoint[
            "model_state_dict"
        ]
    )

    resnet.to(device)


    image_transform = transforms.Compose([
        transforms.Resize(
            (224, 224)
        ),

        transforms.ToTensor(),

        transforms.Normalize(
            mean=[
                0.485,
                0.456,
                0.406
            ],

            std=[
                0.229,
                0.224,
                0.225
            ]
        )
    ])


    # --------------------------------------------------------
    # Export VALIDATION and TEST
    # --------------------------------------------------------

    for split in [
        "validation",
        "test"
    ]:

        print(
            "\n" + "=" * 70
        )

        print(
            split.upper()
        )

        print("=" * 70)

        dataframe = pd.read_parquet(
            DATA_ROOT
            / f"{split}.parquet"
        )

        export_roberta(
            dataframe,
            split,
            roberta,
            tokenizer,
            device
        )

        export_resnet(
            dataframe,
            split,
            resnet,
            image_transform,
            device
        )


    print(
        "\nBaseline probability "
        "export complete."
    )


# END REGISTERED SOURCE BLOCK


In [38]:
%%project_source multimodal-fake-news-detection/scripts/export_baseline_probabilities.py 2
if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


### 5.6 Evaluate late fusion

Join model predictions one-to-one, check labels, search weights using validation macro F1, freeze alpha and evaluate test predictions.

**Source:** `multimodal-fake-news-detection/scripts/evaluate_late_fusion.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `sklearn`  
**Top-level components:** `compute_metrics`, `load_pair`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/baseline_probabilities`
- `results/metrics/late_probability_fusion`

The following cells contain the complete source; Run All registers it for inspection/export.

In [39]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_late_fusion.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd

from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
    confusion_matrix,
)


INPUT_ROOT = Path(
    "results/metrics/baseline_probabilities"
)

OUTPUT_ROOT = Path(
    "results/metrics/late_probability_fusion"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


def compute_metrics(
    labels,
    probabilities
):

    predictions = (
        probabilities >= 0.5
    ).astype(int)

    return {
        "accuracy": float(
            accuracy_score(
                labels,
                predictions
            )
        ),

        "precision": float(
            precision_score(
                labels,
                predictions,
                zero_division=0
            )
        ),

        "recall": float(
            recall_score(
                labels,
                predictions,
                zero_division=0
            )
        ),

        "f1": float(
            f1_score(
                labels,
                predictions,
                zero_division=0
            )
        ),

        "f1_macro": float(
            f1_score(
                labels,
                predictions,
                average="macro",
                zero_division=0
            )
        ),

        "roc_auc": float(
            roc_auc_score(
                labels,
                probabilities
            )
        ),

        "pr_auc": float(
            average_precision_score(
                labels,
                probabilities
            )
        ),

        "confusion_matrix":
            confusion_matrix(
                labels,
                predictions
            ).tolist(),
    }


def load_pair(split):

    roberta = pd.read_csv(
        INPUT_ROOT
        / f"roberta_{split}.csv"
    )

    resnet = pd.read_csv(
        INPUT_ROOT
        / f"resnet_{split}.csv"
    )

    merged = roberta.merge(
        resnet,
        on="id",
        suffixes=(
            "_text",
            "_image"
        ),
        validate="one_to_one"
    )

    if not np.array_equal(
        merged["label_text"],
        merged["label_image"]
    ):

        raise ValueError(
            f"{split}: label mismatch."
        )

    return merged


validation = load_pair(
    "validation"
)

test = load_pair(
    "test"
)


print("=" * 70)
print("LATE PROBABILITY FUSION")
print("=" * 70)

print(
    f"\nValidation samples: "
    f"{len(validation):,}"
)

print(
    f"Test samples:       "
    f"{len(test):,}"
)


# END REGISTERED SOURCE BLOCK


In [40]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_late_fusion.py 1
validation_labels = (
    validation["label_text"]
    .to_numpy()
)

validation_text = (
    validation[
        "probability_class_1_text"
    ]
    .to_numpy()
)

validation_image = (
    validation[
        "probability_class_1_image"
    ]
    .to_numpy()
)


# ------------------------------------------------------------
# Tune alpha ONLY on validation data.
#
# alpha = 1.0 -> text only
# alpha = 0.0 -> image only
# ------------------------------------------------------------

grid_results = []

best_alpha = None
best_macro_f1 = -1.0


for alpha in np.arange(
    0.0,
    1.0001,
    0.05
):

    fused_probability = (
        alpha
        * validation_text
        +
        (1.0 - alpha)
        * validation_image
    )

    metrics = compute_metrics(
        validation_labels,
        fused_probability
    )

    grid_results.append({
        "alpha_text":
            float(round(alpha, 2)),

        "alpha_image":
            float(
                round(
                    1.0 - alpha,
                    2
                )
            ),

        **{
            key: value
            for key, value
            in metrics.items()
            if key !=
            "confusion_matrix"
        }
    })


    current_macro_f1 = (
        metrics["f1_macro"]
    )


    if (
        current_macro_f1
        > best_macro_f1
    ):

        best_macro_f1 = (
            current_macro_f1
        )

        best_alpha = float(
            round(alpha, 2)
        )


grid_df = pd.DataFrame(
    grid_results
)

grid_df.to_csv(
    OUTPUT_ROOT
    / "validation_alpha_search.csv",
    index=False
)


print(
    f"\nBest validation alpha "
    f"(text): {best_alpha:.2f}"
)

print(
    f"Image weight: "
    f"{1.0 - best_alpha:.2f}"
)

print(
    f"Best validation macro F1: "
    f"{best_macro_f1:.4f}"
)


best_validation_probability = (
    best_alpha
    * validation_text
    +
    (1.0 - best_alpha)
    * validation_image
)


validation_metrics = (
    compute_metrics(
        validation_labels,
        best_validation_probability
    )
)


print(
    "\nValidation metrics "
    "at selected alpha:"
)

for key, value in (
    validation_metrics.items()
):

    if key == "confusion_matrix":
        continue

    print(
        f"{key:12s}: "
        f"{value:.4f}"
    )


print(
    "Confusion matrix:"
)

print(
    np.array(
        validation_metrics[
            "confusion_matrix"
        ]
    )
)


# ------------------------------------------------------------
# Freeze alpha.
# Evaluate TEST exactly once.
# ------------------------------------------------------------

# END REGISTERED SOURCE BLOCK


In [41]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_late_fusion.py 2
test_labels = (
    test["label_text"]
    .to_numpy()
)

test_text = (
    test[
        "probability_class_1_text"
    ]
    .to_numpy()
)

test_image = (
    test[
        "probability_class_1_image"
    ]
    .to_numpy()
)


test_probability = (
    best_alpha
    * test_text
    +
    (1.0 - best_alpha)
    * test_image
)


test_metrics = compute_metrics(
    test_labels,
    test_probability
)


print("\n" + "=" * 70)
print("TEST RESULTS")
print("=" * 70)


for key, value in (
    test_metrics.items()
):

    if key == "confusion_matrix":
        continue

    print(
        f"{key:12s}: "
        f"{value:.4f}"
    )


print(
    "\nConfusion matrix:"
)

print(
    np.array(
        test_metrics[
            "confusion_matrix"
        ]
    )
)


test_predictions = (
    test_probability >= 0.5
).astype(int)


pd.DataFrame({
    "id":
        test["id"],

    "label":
        test_labels,

    "probability_text":
        test_text,

    "probability_image":
        test_image,

    "probability_fused":
        test_probability,

    "prediction":
        test_predictions,
}).to_csv(
    OUTPUT_ROOT
    / "test_predictions.csv",
    index=False
)


with (
    OUTPUT_ROOT
    / "results.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        {
            "selected_alpha_text":
                best_alpha,

            "selected_alpha_image":
                1.0 - best_alpha,

            "selection_metric":
                "validation_macro_f1",

            "validation":
                validation_metrics,

            "test":
                test_metrics,
        },

        f,
        indent=2
    )


print(
    "\nResults saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


<a id="diagnostics"></a>
## 6. Development diagnostics and explainability

These original diagnostic scripts consume development artifacts. Final-holdout statistics are also produced separately in the next section.

### 6.1 Compare fusion vs roberta

Compare paired development predictions using the implemented statistical tests and bootstrap calculations.

**Source:** `multimodal-fake-news-detection/scripts/compare_fusion_vs_roberta.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `scipy`, `sklearn`  
**Top-level components:** `calculate_metrics`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/baseline_probabilities`
- `results/metrics/late_probability_fusion`
- `results/metrics/statistical_comparison`

The following cells contain the complete source; Run All registers it for inspection/export.

In [42]:
%%project_source multimodal-fake-news-detection/scripts/compare_fusion_vs_roberta.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd

from scipy.stats import binomtest

from sklearn.metrics import (
    accuracy_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
)


SEED = 42
N_BOOTSTRAPS = 5000

BASELINE_ROOT = Path(
    "results/metrics/baseline_probabilities"
)

FUSION_ROOT = Path(
    "results/metrics/late_probability_fusion"
)

OUTPUT_ROOT = Path(
    "results/metrics/statistical_comparison"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


# ============================================================
# Load paired predictions
# ============================================================

roberta = pd.read_csv(
    BASELINE_ROOT / "roberta_test.csv"
)

fusion = pd.read_csv(
    FUSION_ROOT / "test_predictions.csv"
)


df = roberta.merge(
    fusion,
    on="id",
    suffixes=("_roberta", "_fusion"),
    validate="one_to_one"
)


if not np.array_equal(
    df["label_roberta"],
    df["label_fusion"]
):
    raise ValueError(
        "Label mismatch between prediction files."
    )


y = df["label_roberta"].to_numpy()

pred_roberta = (
    df["prediction_roberta"]
    .to_numpy()
)

pred_fusion = (
    df["prediction_fusion"]
    .to_numpy()
)

prob_roberta = (
    df["probability_class_1"]
    .to_numpy()
)

prob_fusion = (
    df["probability_fused"]
    .to_numpy()
)


print("=" * 70)
print("LATE FUSION VS ROBERTA")
print("=" * 70)

print(f"\nPaired test samples: {len(df):,}")


# ============================================================
# McNemar exact test
# ============================================================

correct_roberta = (
    pred_roberta == y
)

correct_fusion = (
    pred_fusion == y
)


# RoBERTa correct, fusion wrong
b = int(
    np.sum(
        correct_roberta
        & ~correct_fusion
    )
)

# RoBERTa wrong, fusion correct
c = int(
    np.sum(
        ~correct_roberta
        & correct_fusion
    )
)


discordant = b + c


if discordant > 0:

    mcnemar = binomtest(
        min(b, c),
        n=discordant,
        p=0.5,
        alternative="two-sided"
    )

    mcnemar_p = float(
        mcnemar.pvalue
    )

else:
    mcnemar_p = 1.0


print("\nMcNemar paired comparison:")
print(
    "RoBERTa correct / Fusion wrong:",
    b
)

print(
    "RoBERTa wrong / Fusion correct:",
    c
)

print(
    "Discordant predictions:",
    discordant
)

# END REGISTERED SOURCE BLOCK


In [43]:
%%project_source multimodal-fake-news-detection/scripts/compare_fusion_vs_roberta.py 1
print(
    f"Exact p-value: {mcnemar_p:.6f}"
)


# ============================================================
# Metric helper
# ============================================================

def calculate_metrics(
    labels,
    predictions,
    probabilities
):

    return {
        "accuracy":
            accuracy_score(
                labels,
                predictions
            ),

        "f1":
            f1_score(
                labels,
                predictions
            ),

        "f1_macro":
            f1_score(
                labels,
                predictions,
                average="macro"
            ),

        "roc_auc":
            roc_auc_score(
                labels,
                probabilities
            ),

        "pr_auc":
            average_precision_score(
                labels,
                probabilities
            ),
    }


roberta_metrics = calculate_metrics(
    y,
    pred_roberta,
    prob_roberta
)

fusion_metrics = calculate_metrics(
    y,
    pred_fusion,
    prob_fusion
)


print("\nObserved metric differences:")
print("(Fusion - RoBERTa)")

for metric in roberta_metrics:

    delta = (
        fusion_metrics[metric]
        - roberta_metrics[metric]
    )

    print(
        f"{metric:12s}: "
        f"{delta:+.4f}"
    )


# ============================================================
# Paired bootstrap
# ============================================================

rng = np.random.default_rng(
    SEED
)

n = len(df)

bootstrap_differences = {
    metric: []
    for metric in roberta_metrics
}


print(
    f"\nRunning {N_BOOTSTRAPS:,} "
    "paired bootstrap samples..."
)


for i in range(N_BOOTSTRAPS):

    indices = rng.integers(
        0,
        n,
        size=n
    )

    y_sample = y[indices]

    # ROC/PR require both labels to appear.
    if len(np.unique(y_sample)) < 2:
        continue

    roberta_sample = (
        calculate_metrics(
            y_sample,
            pred_roberta[indices],
            prob_roberta[indices]
        )
    )

    fusion_sample = (
        calculate_metrics(
            y_sample,
            pred_fusion[indices],
            prob_fusion[indices]
        )
    )

    for metric in (
        bootstrap_differences
    ):

        bootstrap_differences[
            metric
        ].append(
            fusion_sample[metric]
            - roberta_sample[metric]
        )


# ============================================================
# Confidence intervals
# ============================================================

confidence_intervals = {}


print("\n95% bootstrap confidence intervals:")
print("(Fusion - RoBERTa)")


for metric, differences in (
    bootstrap_differences.items()
):

    values = np.asarray(
        differences
    )

    lower = float(
        np.percentile(
            values,
            2.5
        )
    )

    upper = float(
        np.percentile(
            values,
            97.5
        )
    )

    observed = float(
        fusion_metrics[metric]
        - roberta_metrics[metric]
    )

    confidence_intervals[
        metric
    ] = {
        "observed_difference":
            observed,

        "ci_95_lower":
            lower,

        "ci_95_upper":
            upper,
    }

    print(
        f"{metric:12s}: "
        f"{observed:+.4f} "
        f"[{lower:+.4f}, {upper:+.4f}]"
    )


# ============================================================
# Save results
# ============================================================

# END REGISTERED SOURCE BLOCK


In [44]:
%%project_source multimodal-fake-news-detection/scripts/compare_fusion_vs_roberta.py 2
results = {
    "comparison":
        "late_probability_fusion_vs_roberta",

    "test_samples":
        int(n),

    "mcnemar": {
        "roberta_correct_fusion_wrong":
            b,

        "roberta_wrong_fusion_correct":
            c,

        "discordant":
            discordant,

        "exact_p_value":
            mcnemar_p,
    },

    "roberta_metrics": {
        key: float(value)
        for key, value
        in roberta_metrics.items()
    },

    "fusion_metrics": {
        key: float(value)
        for key, value
        in fusion_metrics.items()
    },

    "bootstrap_samples":
        N_BOOTSTRAPS,

    "confidence_intervals":
        confidence_intervals,
}


with (
    OUTPUT_ROOT / "results.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        results,
        f,
        indent=2
    )


print(
    "\nResults saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


### 6.2 Analyse calibration

Measure whether predictive probabilities agree with empirical outcomes, using Brier score, log loss and calibration summaries.

**Source:** `multimodal-fake-news-detection/scripts/analyse_calibration.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `sklearn`  
**Top-level components:** `expected_calibration_error`, `model_calibration`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/baseline_probabilities`
- `results/metrics/late_probability_fusion`
- `results/metrics/calibration_analysis`

The following cells contain the complete source; Run All registers it for inspection/export.

In [45]:
%%project_source multimodal-fake-news-detection/scripts/analyse_calibration.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd

from sklearn.metrics import (
    brier_score_loss,
    log_loss,
)


PROB_ROOT = Path(
    "results/metrics/baseline_probabilities"
)

FUSION_ROOT = Path(
    "results/metrics/late_probability_fusion"
)

OUTPUT_ROOT = Path(
    "results/metrics/calibration_analysis"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


N_BINS = 10


def expected_calibration_error(
    labels,
    probabilities,
    n_bins=10
):

    probabilities = np.asarray(
        probabilities
    )

    labels = np.asarray(
        labels
    )

    predictions = (
        probabilities >= 0.5
    ).astype(int)

    confidence = np.maximum(
        probabilities,
        1.0 - probabilities
    )

    correctness = (
        predictions == labels
    ).astype(float)

    bin_edges = np.linspace(
        0.5,
        1.0,
        n_bins + 1
    )

    ece = 0.0
    rows = []

    for i in range(n_bins):

        lower = bin_edges[i]
        upper = bin_edges[i + 1]

        if i == n_bins - 1:
            mask = (
                (confidence >= lower)
                & (confidence <= upper)
            )
        else:
            mask = (
                (confidence >= lower)
                & (confidence < upper)
            )

        count = int(mask.sum())

        if count == 0:
            rows.append({
                "bin_lower": lower,
                "bin_upper": upper,
                "count": 0,
                "mean_confidence": None,
                "accuracy": None,
                "gap": None,
            })

            continue

        mean_confidence = float(
            confidence[mask].mean()
        )

        accuracy = float(
            correctness[mask].mean()
        )

        gap = abs(
            accuracy - mean_confidence
        )

        ece += (
            count / len(labels)
        ) * gap

        rows.append({
            "bin_lower": float(lower),
            "bin_upper": float(upper),
            "count": count,
            "mean_confidence":
                mean_confidence,
            "accuracy":
                accuracy,
            "gap":
                float(gap),
        })

    return float(ece), rows


def model_calibration(
    name,
    labels,
    probabilities
):

    probabilities = np.clip(
        np.asarray(probabilities),
        1e-7,
        1 - 1e-7
    )

    ece, bins = (
        expected_calibration_error(
            labels,
            probabilities,
            N_BINS
        )
    )

    result = {
        "model": name,

        "brier_score":
            float(
                brier_score_loss(
                    labels,
                    probabilities
                )
            ),

        "log_loss":
            float(
                log_loss(
                    labels,
                    probabilities
                )
            ),

        "ece":
            ece,

        "mean_probability_class_1":
            float(
                probabilities.mean()
            ),

        "mean_confidence":
            float(
                np.maximum(
                    probabilities,
                    1 - probabilities
                ).mean()
            ),
    }

    return result, bins


# END REGISTERED SOURCE BLOCK


In [46]:
%%project_source multimodal-fake-news-detection/scripts/analyse_calibration.py 1
roberta = pd.read_csv(
    PROB_ROOT / "roberta_test.csv"
)

resnet = pd.read_csv(
    PROB_ROOT / "resnet_test.csv"
)

fusion = pd.read_csv(
    FUSION_ROOT / "test_predictions.csv"
)


df = (
    roberta[
        [
            "id",
            "label",
            "probability_class_1"
        ]
    ]
    .rename(
        columns={
            "probability_class_1":
                "probability_roberta"
        }
    )
    .merge(
        resnet[
            [
                "id",
                "probability_class_1"
            ]
        ].rename(
            columns={
                "probability_class_1":
                    "probability_resnet"
            }
        ),
        on="id",
        validate="one_to_one"
    )
    .merge(
        fusion[
            [
                "id",
                "probability_fused"
            ]
        ],
        on="id",
        validate="one_to_one"
    )
)


labels = (
    df["label"]
    .to_numpy()
)


models = {
    "roberta":
        df[
            "probability_roberta"
        ].to_numpy(),

    "resnet":
        df[
            "probability_resnet"
        ].to_numpy(),

    "late_fusion":
        df[
            "probability_fused"
        ].to_numpy(),
}


summary = []
all_bins = {}


print("=" * 70)
print("MODEL CALIBRATION ANALYSIS")
print("=" * 70)

print(
    f"\nTest samples: {len(df):,}"
)


for name, probabilities in (
    models.items()
):

    result, bins = (
        model_calibration(
            name,
            labels,
            probabilities
        )
    )

    summary.append(
        result
    )

    all_bins[name] = bins

    print(
        "\n" + name.upper()
    )

    print(
        "-" * len(name)
    )

    print(
        f"Brier score : "
        f"{result['brier_score']:.4f}"
    )

    print(
        f"Log loss    : "
        f"{result['log_loss']:.4f}"
    )

    print(
        f"ECE         : "
        f"{result['ece']:.4f}"
    )

    print(
        f"Mean conf.  : "
        f"{result['mean_confidence']:.4f}"
    )


summary_df = pd.DataFrame(
    summary
)

summary_df.to_csv(
    OUTPUT_ROOT
    / "calibration_summary.csv",
    index=False
)


for model, bins in (
    all_bins.items()
):

    pd.DataFrame(
        bins
    ).to_csv(
        OUTPUT_ROOT
        / f"{model}_calibration_bins.csv",
        index=False
    )


# END REGISTERED SOURCE BLOCK


In [47]:
%%project_source multimodal-fake-news-detection/scripts/analyse_calibration.py 2
with (
    OUTPUT_ROOT
    / "results.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        {
            "n_bins":
                N_BINS,

            "test_samples":
                int(len(df)),

            "models":
                summary,
        },
        f,
        indent=2
    )


print(
    "\n" + "=" * 70
)

print(
    "SUMMARY"
)

print("=" * 70)

print(
    summary_df[
        [
            "model",
            "brier_score",
            "log_loss",
            "ece",
            "mean_confidence",
        ]
    ].to_string(
        index=False,
        float_format=lambda x:
            f"{x:.4f}"
    )
)

print(
    "\nLower Brier, log loss, "
    "and ECE indicate better calibration."
)

print(
    "\nResults saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


### 6.3 Analyse missing modality

Study the implemented missing-modality conditions and fallback behaviour; distinguish simulated removal from naturally absent images.

**Source:** `multimodal-fake-news-detection/scripts/analyse_missing_modality.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `sklearn`  
**Top-level components:** `metrics`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/baseline_probabilities`
- `results/metrics/missing_modality_robustness`

The following cells contain the complete source; Run All registers it for inspection/export.

In [48]:
%%project_source multimodal-fake-news-detection/scripts/analyse_missing_modality.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd

from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
)


INPUT_ROOT = Path(
    "results/metrics/baseline_probabilities"
)

OUTPUT_ROOT = Path(
    "results/metrics/missing_modality_robustness"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


ALPHA_TEXT = 0.45
ALPHA_IMAGE = 0.55

THRESHOLD = 0.5


def metrics(
    labels,
    probabilities
):

    predictions = (
        probabilities >= THRESHOLD
    ).astype(int)

    return {
        "accuracy":
            float(
                accuracy_score(
                    labels,
                    predictions
                )
            ),

        "precision":
            float(
                precision_score(
                    labels,
                    predictions,
                    zero_division=0
                )
            ),

        "recall":
            float(
                recall_score(
                    labels,
                    predictions,
                    zero_division=0
                )
            ),

        "f1":
            float(
                f1_score(
                    labels,
                    predictions,
                    zero_division=0
                )
            ),

        "f1_macro":
            float(
                f1_score(
                    labels,
                    predictions,
                    average="macro",
                    zero_division=0
                )
            ),

        "roc_auc":
            float(
                roc_auc_score(
                    labels,
                    probabilities
                )
            ),

        "pr_auc":
            float(
                average_precision_score(
                    labels,
                    probabilities
                )
            ),
    }


# ============================================================
# VALIDATION ONLY
# ============================================================

text = pd.read_csv(
    INPUT_ROOT
    / "roberta_validation.csv"
)

image = pd.read_csv(
    INPUT_ROOT
    / "resnet_validation.csv"
)


df = text.merge(
    image,
    on="id",
    suffixes=(
        "_text",
        "_image"
    ),
    validate="one_to_one"
)


if not np.array_equal(
    df["label_text"],
    df["label_image"]
):

    raise ValueError(
        "Validation labels do not match."
    )


labels = (
    df["label_text"]
    .to_numpy()
)

p_text = (
    df[
        "probability_class_1_text"
    ]
    .to_numpy()
)

p_image = (
    df[
        "probability_class_1_image"
    ]
    .to_numpy()
)


# ============================================================
# Scenarios
# ============================================================

# END REGISTERED SOURCE BLOCK


In [49]:
%%project_source multimodal-fake-news-detection/scripts/analyse_missing_modality.py 1
scenarios = {}


# Full multimodal model
scenarios["normal_late_fusion"] = (
    ALPHA_TEXT
    * p_text
    +
    ALPHA_IMAGE
    * p_image
)


# Explicit fallback strategies
scenarios["missing_image_text_fallback"] = (
    p_text
)

scenarios["missing_text_image_fallback"] = (
    p_image
)


# Naive neutral-imputation strategies
scenarios["missing_image_neutral"] = (
    ALPHA_TEXT
    * p_text
    +
    ALPHA_IMAGE
    * 0.5
)

scenarios["missing_text_neutral"] = (
    ALPHA_TEXT
    * 0.5
    +
    ALPHA_IMAGE
    * p_image
)


# ============================================================
# Evaluate
# ============================================================

results = []


print("=" * 70)
print("MISSING-MODALITY ROBUSTNESS")
print("=" * 70)

print(
    f"\nValidation samples: "
    f"{len(df):,}"
)

print(
    "\nTEST SET IS NOT USED."
)


for name, probability in (
    scenarios.items()
):

    result = metrics(
        labels,
        probability
    )

    result["scenario"] = name

    results.append(
        result
    )


    print(
        "\n" + name.upper()
    )

    print(
        "-" * len(name)
    )

    for metric, value in (
        result.items()
    ):

        if metric == "scenario":
            continue

        print(
            f"{metric:12s}: "
            f"{value:.4f}"
        )


results_df = pd.DataFrame(
    results
)


baseline_macro = float(
    results_df.loc[
        results_df["scenario"]
        == "normal_late_fusion",
        "f1_macro"
    ].iloc[0]
)


results_df[
    "macro_f1_change_vs_full"
] = (
    results_df["f1_macro"]
    - baseline_macro
)


results_df.to_csv(
    OUTPUT_ROOT
    / "robustness_results.csv",
    index=False
)


with (
    OUTPUT_ROOT
    / "results.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        {
            "dataset_split":
                "validation",

            "test_used":
                False,

            "alpha_text":
                ALPHA_TEXT,

            "alpha_image":
                ALPHA_IMAGE,

            "results":
                results_df
                .to_dict(
                    orient="records"
                ),
        },
        f,
        indent=2
    )


# END REGISTERED SOURCE BLOCK


In [50]:
%%project_source multimodal-fake-news-detection/scripts/analyse_missing_modality.py 2
print(
    "\n" + "=" * 70
)

print(
    "SUMMARY"
)

print("=" * 70)

print(
    results_df[
        [
            "scenario",
            "accuracy",
            "f1_macro",
            "roc_auc",
            "pr_auc",
            "macro_f1_change_vs_full",
        ]
    ].to_string(
        index=False,
        float_format=lambda x:
            f"{x:.4f}"
    )
)


print(
    "\nResults saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


### 6.4 Analyse model errors

Identify agreement/disagreement patterns and examples where one modality helps or hurts.

**Source:** `multimodal-fake-news-detection/scripts/analyse_model_errors.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/baseline_probabilities`
- `results/metrics/late_probability_fusion`
- `data/processed/fakeddit/development_clean/test.parquet`
- `results/metrics/error_analysis`

The following cells contain the complete source; Run All registers it for inspection/export.

In [51]:
%%project_source multimodal-fake-news-detection/scripts/analyse_model_errors.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd


PROB_ROOT = Path(
    "results/metrics/baseline_probabilities"
)

FUSION_ROOT = Path(
    "results/metrics/late_probability_fusion"
)

DATA_PATH = Path(
    "data/processed/fakeddit/development_clean/test.parquet"
)

OUTPUT_ROOT = Path(
    "results/metrics/error_analysis"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


roberta = pd.read_csv(
    PROB_ROOT / "roberta_test.csv"
)

resnet = pd.read_csv(
    PROB_ROOT / "resnet_test.csv"
)

fusion = pd.read_csv(
    FUSION_ROOT / "test_predictions.csv"
)

data = pd.read_parquet(
    DATA_PATH
)


# ------------------------------------------------------------
# Standardise IDs
# ------------------------------------------------------------

for frame in [
    roberta,
    resnet,
    fusion,
    data
]:
    frame["id"] = (
        frame["id"]
        .astype(str)
    )


# ------------------------------------------------------------
# Rename model outputs
# ------------------------------------------------------------

roberta = roberta.rename(
    columns={
        "prediction":
            "prediction_roberta",

        "probability_class_1":
            "probability_roberta",
    }
)

resnet = resnet.rename(
    columns={
        "prediction":
            "prediction_resnet",

        "probability_class_1":
            "probability_resnet",
    }
)

fusion = fusion.rename(
    columns={
        "prediction":
            "prediction_fusion",
    }
)


# ------------------------------------------------------------
# Merge paired results
# ------------------------------------------------------------

df = (
    data
    .merge(
        roberta[
            [
                "id",
                "prediction_roberta",
                "probability_roberta",
            ]
        ],
        on="id",
        validate="one_to_one"
    )
    .merge(
        resnet[
            [
                "id",
                "prediction_resnet",
                "probability_resnet",
            ]
        ],
        on="id",
        validate="one_to_one"
    )
    .merge(
        fusion[
            [
                "id",
                "prediction_fusion",
                "probability_fused",
            ]
        ],
        on="id",
        validate="one_to_one"
    )
)


df["roberta_correct"] = (
    df["prediction_roberta"]
    == df["label"]
)

df["resnet_correct"] = (
    df["prediction_resnet"]
    == df["label"]
)

df["fusion_correct"] = (
    df["prediction_fusion"]
    == df["label"]
)


# ------------------------------------------------------------
# Pairwise categories
# ------------------------------------------------------------

conditions = [
    (
        df["roberta_correct"]
        & df["fusion_correct"]
    ),

    (
        ~df["roberta_correct"]
        & df["fusion_correct"]
    ),

    (
        df["roberta_correct"]
        & ~df["fusion_correct"]
    ),

    (
        ~df["roberta_correct"]
        & ~df["fusion_correct"]
    ),
]

# END REGISTERED SOURCE BLOCK


In [52]:
%%project_source multimodal-fake-news-detection/scripts/analyse_model_errors.py 1
categories = [
    "both_correct",
    "fusion_only_correct",
    "roberta_only_correct",
    "both_wrong",
]

df["comparison_group"] = np.select(
    conditions,
    categories,
    default="unknown"
)


# ------------------------------------------------------------
# Basic counts
# ------------------------------------------------------------

counts = (
    df["comparison_group"]
    .value_counts()
    .to_dict()
)

print("=" * 70)
print("ERROR / COMPLEMENTARITY ANALYSIS")
print("=" * 70)

print("\nRoBERTa vs Fusion groups:")

for group in categories:
    print(
        f"{group:22s}: "
        f"{counts.get(group, 0):,}"
    )


# ------------------------------------------------------------
# Recovered cases
# ------------------------------------------------------------

recovered = df[
    df["comparison_group"]
    == "fusion_only_correct"
].copy()

lost = df[
    df["comparison_group"]
    == "roberta_only_correct"
].copy()


print("\nFusion recovered cases:")
print(
    f"Total: {len(recovered):,}"
)

print("\nRecovered cases by true label:")
print(
    recovered["label"]
    .value_counts()
    .sort_index()
)


resnet_correct_recovered = int(
    recovered[
        "resnet_correct"
    ].sum()
)


print(
    "\nAmong recovered cases, "
    "ResNet was independently correct:"
)

print(
    f"{resnet_correct_recovered:,} "
    f"/ {len(recovered):,} "
    f"("
    f"{resnet_correct_recovered / len(recovered):.1%}"
    f")"
)


print("\nFusion-lost cases:")
print(
    f"Total: {len(lost):,}"
)

print("\nLost cases by true label:")
print(
    lost["label"]
    .value_counts()
    .sort_index()
)


# ------------------------------------------------------------
# Model agreement
# ------------------------------------------------------------

agreement = (
    df["prediction_roberta"]
    == df["prediction_resnet"]
)

print(
    "\nRoBERTa / ResNet prediction agreement:"
)

print(
    f"{agreement.mean():.1%}"
)


disagreement = df[
    ~agreement
].copy()

print(
    "Samples where modalities disagree:",
    len(disagreement)
)

print(
    "\nWhen RoBERTa and ResNet disagree:"
)

print(
    "RoBERTa correct:",
    int(
        disagreement[
            "roberta_correct"
        ].sum()
    )
)

print(
    "ResNet correct:",
    int(
        disagreement[
            "resnet_correct"
        ].sum()
    )
)

print(
    "Fusion correct:",
    int(
        disagreement[
            "fusion_correct"
        ].sum()
    )
)


# ------------------------------------------------------------
# Text length
# ------------------------------------------------------------

# END REGISTERED SOURCE BLOCK


In [53]:
%%project_source multimodal-fake-news-detection/scripts/analyse_model_errors.py 2
if "text_length_words" in df.columns:
    text_length = "text_length_words"
else:
    df["derived_text_words"] = (
        df["text"]
        .fillna("")
        .astype(str)
        .str.split()
        .str.len()
    )

    text_length = (
        "derived_text_words"
    )


print("\nMean text length by group:")

print(
    df.groupby(
        "comparison_group"
    )[text_length]
    .mean()
    .reindex(categories)
)


# ------------------------------------------------------------
# Probability shifts
# ------------------------------------------------------------

df[
    "fusion_minus_roberta_probability"
] = (
    df["probability_fused"]
    - df["probability_roberta"]
)


print(
    "\nMean probability shift "
    "(Fusion - RoBERTa) by group:"
)

print(
    df.groupby(
        "comparison_group"
    )[
        "fusion_minus_roberta_probability"
    ]
    .mean()
    .reindex(categories)
)


# ------------------------------------------------------------
# Save detailed data
# ------------------------------------------------------------

df.to_csv(
    OUTPUT_ROOT
    / "paired_test_error_analysis.csv",
    index=False
)

recovered.to_csv(
    OUTPUT_ROOT
    / "fusion_recovered_cases.csv",
    index=False
)

lost.to_csv(
    OUTPUT_ROOT
    / "fusion_lost_cases.csv",
    index=False
)


summary = {
    "test_samples":
        int(len(df)),

    "groups": {
        key: int(value)
        for key, value
        in counts.items()
    },

    "fusion_recovered":
        int(len(recovered)),

    "fusion_lost":
        int(len(lost)),

    "resnet_correct_among_recovered":
        resnet_correct_recovered,

    "resnet_correct_among_recovered_rate":
        float(
            resnet_correct_recovered
            / len(recovered)
        ),

    "roberta_resnet_agreement":
        float(
            agreement.mean()
        ),

    "modality_disagreement_samples":
        int(len(disagreement)),

    "when_modalities_disagree": {
        "roberta_correct":
            int(
                disagreement[
                    "roberta_correct"
                ].sum()
            ),

        "resnet_correct":
            int(
                disagreement[
                    "resnet_correct"
                ].sum()
            ),

        "fusion_correct":
            int(
                disagreement[
                    "fusion_correct"
                ].sum()
            ),
    },
}


with (
    OUTPUT_ROOT / "summary.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        summary,
        f,
        indent=2
    )


print(
    "\nResults saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


### 6.5 Generate roberta shap cases

Generate selected text attributions from the saved model. These are explanations of model behaviour, not proof of factual validity.

**Source:** `multimodal-fake-news-detection/scripts/generate_roberta_shap_cases.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`, `shap`, `torch`, `transformers`  
**Top-level components:** `predict_proba`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `checkpoints/roberta_baseline`
- `results/gradcam/gradcam_case_summary.csv`
- `results/shap`

The following cells contain the complete source; Run All registers it for inspection/export.

In [54]:
%%project_source multimodal-fake-news-detection/scripts/generate_roberta_shap_cases.py 0
from pathlib import Path
import json

import numpy as np
import pandas as pd
import torch
import shap

from transformers import (
    AutoTokenizer,
    AutoModelForSequenceClassification,
)


CHECKPOINT_PATH = Path(
    "checkpoints/roberta_baseline"
)

CASE_PATH = Path(
    "results/gradcam/gradcam_case_summary.csv"
)

OUTPUT_ROOT = Path(
    "results/shap"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


MAX_LENGTH = 64
MAX_EVALS = 128
BATCH_SIZE = 32


device = torch.device(
    "cuda"
    if torch.cuda.is_available()
    else "cpu"
)


print("=" * 70)
print("ROBERTA SHAP TEXT ATTRIBUTION")
print("=" * 70)

print(
    f"\nDevice: {device}"
)

if device.type == "cuda":

    print(
        "GPU:",
        torch.cuda.get_device_name(0)
    )


# ============================================================
# Load fine-tuned RoBERTa
# ============================================================

print(
    "\nLoading RoBERTa checkpoint..."
)

tokenizer = (
    AutoTokenizer
    .from_pretrained(
        CHECKPOINT_PATH
    )
)

model = (
    AutoModelForSequenceClassification
    .from_pretrained(
        CHECKPOINT_PATH
    )
)

model.to(device)
model.eval()


# ============================================================
# Prediction function used by SHAP
# ============================================================

def predict_proba(texts):

    texts = [
        str(text)
        for text in texts
    ]

    encoded = tokenizer(
        texts,
        padding=True,
        truncation=True,
        max_length=MAX_LENGTH,
        return_tensors="pt"
    )

    encoded = {
        key: value.to(device)
        for key, value
        in encoded.items()
    }

    with torch.no_grad():

        logits = model(
            **encoded
        ).logits

        probabilities = torch.softmax(
            logits,
            dim=1
        )

    return (
        probabilities
        .cpu()
        .numpy()
    )


# ============================================================
# SHAP explainer
# ============================================================

masker = shap.maskers.Text(
    tokenizer
)

explainer = shap.Explainer(
    predict_proba,
    masker,
    algorithm="partition",
    output_names=[
        "class_0",
        "class_1",
    ]
)


# ============================================================
# Load same 32 cases as Grad-CAM
# ============================================================

cases = pd.read_csv(
    CASE_PATH
)

print(
    f"\nCases: {len(cases):,}"
)


# END REGISTERED SOURCE BLOCK


In [55]:
%%project_source multimodal-fake-news-detection/scripts/generate_roberta_shap_cases.py 1
all_token_rows = []
case_summaries = []


for index, row in cases.iterrows():

    sample_id = str(
        row["id"]
    )

    text = str(
        row["text"]
    )

    expected_prediction = int(
        row["prediction_roberta"]
    )


    print(
        "\n" + "=" * 70
    )

    print(
        f"{index + 1}/{len(cases)} "
        f"{sample_id}"
    )

    print(
        f"Group: "
        f"{row['comparison_group']}"
    )

    print(
        f"Text: {text}"
    )


    # --------------------------------------------------------
    # Verify current model prediction
    # --------------------------------------------------------

    probability = predict_proba(
        [text]
    )[0]

    predicted_class = int(
        np.argmax(
            probability
        )
    )


    print(
        "Probability class 0:",
        f"{probability[0]:.4f}"
    )

    print(
        "Probability class 1:",
        f"{probability[1]:.4f}"
    )

    print(
        "Predicted class:",
        predicted_class
    )


    if (
        predicted_class
        != expected_prediction
    ):

        print(
            "WARNING: prediction differs "
            "from stored evaluation output."
        )


    # --------------------------------------------------------
    # SHAP explanation
    #
    # We explain the class actually predicted
    # by RoBERTa.
    # --------------------------------------------------------

    explanation = explainer(
        [text],
        max_evals=MAX_EVALS,
        batch_size=BATCH_SIZE
    )


    tokens = list(
        explanation.data[0]
    )

    values = (
        explanation.values[
            0,
            :,
            predicted_class
        ]
    )


    # --------------------------------------------------------
    # Save token attributions
    # --------------------------------------------------------

    token_rows = []


    for token, value in zip(
        tokens,
        values
    ):

        cleaned_token = str(
            token
        )

        attribution = float(
            value
        )


        token_row = {
            "id":
                sample_id,

            "comparison_group":
                row[
                    "comparison_group"
                ],

            "label":
                int(
                    row["label"]
                ),

            "predicted_class":
                predicted_class,

            "token":
                cleaned_token,

            "shap_value":
                attribution,

            "absolute_shap":
                abs(attribution),
        }


        token_rows.append(
            token_row
        )

        all_token_rows.append(
            token_row
        )


    token_df = pd.DataFrame(
        token_rows
    )


    token_df.to_csv(
        OUTPUT_ROOT
        / f"{sample_id}_tokens.csv",
        index=False
    )


    # --------------------------------------------------------
    # Top supportive/opposing tokens
    # --------------------------------------------------------

    meaningful = token_df[
        token_df["token"]
        .astype(str)
        .str.strip()
        .ne("")
    ].copy()


    supportive = (
        meaningful
        .sort_values(
            "shap_value",
            ascending=False
        )
        .head(5)
    )


    opposing = (
        meaningful
        .sort_values(
            "shap_value",
            ascending=True
        )
        .head(5)
    )


    supportive_text = [
        {
            "token":
                str(r["token"]),

            "value":
                float(
                    r["shap_value"]
                ),
        }

        for _, r
        in supportive.iterrows()
    ]


    opposing_text = [
        {
            "token":
                str(r["token"]),

            "value":
                float(
                    r["shap_value"]
                ),
        }

        for _, r
        in opposing.iterrows()
    ]


    print(
        "\nTop tokens supporting "
        f"class {predicted_class}:"
    )

    for item in supportive_text:

        print(
            f"  {item['token']!r}: "
            f"{item['value']:+.4f}"
        )


    print(
        "\nTop tokens opposing "
        f"class {predicted_class}:"
    )

    for item in opposing_text:

        print(
            f"  {item['token']!r}: "
            f"{item['value']:+.4f}"
        )


    case_summaries.append({
        "id":
            sample_id,

        "comparison_group":
            row[
                "comparison_group"
            ],

        "text":
            text,

        "label":
            int(
                row["label"]
            ),

        "prediction_roberta":
            expected_prediction,

        "shap_predicted_class":
            predicted_class,

        "probability_class_0":
            float(
                probability[0]
            ),

        "probability_class_1":
            float(
                probability[1]
            ),

        "top_supportive_tokens":
            json.dumps(
                supportive_text
            ),

        "top_opposing_tokens":
            json.dumps(
                opposing_text
            ),
    })


# ============================================================
# Save consolidated outputs
# ============================================================

# END REGISTERED SOURCE BLOCK


In [56]:
%%project_source multimodal-fake-news-detection/scripts/generate_roberta_shap_cases.py 2
pd.DataFrame(
    all_token_rows
).to_csv(
    OUTPUT_ROOT
    / "all_token_attributions.csv",
    index=False
)


pd.DataFrame(
    case_summaries
).to_csv(
    OUTPUT_ROOT
    / "shap_case_summary.csv",
    index=False
)


with (
    OUTPUT_ROOT
    / "metadata.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        {
            "method":
                "SHAP Partition Explainer",

            "model":
                "fine-tuned roberta-base",

            "cases":
                int(len(cases)),

            "max_length":
                MAX_LENGTH,

            "max_evals":
                MAX_EVALS,

            "explained_output":
                "RoBERTa predicted class",

            "interpretation":
                (
                    "Positive SHAP values support "
                    "the predicted class; negative "
                    "values oppose the predicted class."
                ),
        },
        f,
        indent=2
    )


print(
    "\n" + "=" * 70
)

print(
    "ROBERTA SHAP COMPLETE"
)

print("=" * 70)

print(
    f"\nExplained {len(cases):,} cases."
)

print(
    "Saved to:",
    OUTPUT_ROOT
)


if __name__ == "__main__":
    pass
# END REGISTERED SOURCE BLOCK


### 6.6 Generate gradcam cases

Generate selected visual activation explanations using the saved image model.

**Source:** `multimodal-fake-news-detection/scripts/generate_gradcam_cases.py`  
**Imported modules:** `PIL`, `numpy`, `pandas`, `pathlib`, `pytorch_grad_cam`, `random`, `torch`, `torchvision`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/metrics/error_analysis/paired_test_error_analysis.csv`
- `checkpoints/resnet50_baseline/best_model.pt`
- `results/gradcam`

The following cells contain the complete source; Run All registers it for inspection/export.

In [57]:
%%project_source multimodal-fake-news-detection/scripts/generate_gradcam_cases.py 0
from pathlib import Path
import random

import numpy as np
import pandas as pd
from PIL import Image
from pytorch_grad_cam.utils.model_targets import (
    ClassifierOutputTarget,
)

import torch
import torch.nn as nn

from torchvision.models import resnet50
from torchvision import transforms

from pytorch_grad_cam import GradCAM
from pytorch_grad_cam.utils.image import (
    show_cam_on_image,
)


SEED = 42
N_PER_GROUP = 8

ERROR_PATH = Path(
    "results/metrics/error_analysis/"
    "paired_test_error_analysis.csv"
)

CHECKPOINT_PATH = Path(
    "checkpoints/resnet50_baseline/best_model.pt"
)

OUTPUT_ROOT = Path(
    "results/gradcam"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


random.seed(SEED)
np.random.seed(SEED)
torch.manual_seed(SEED)


device = torch.device(
    "cuda"
    if torch.cuda.is_available()
    else "cpu"
)


# ============================================================
# Load ResNet
# ============================================================

model = resnet50(
    weights=None
)

features = model.fc.in_features

model.fc = nn.Linear(
    features,
    2
)


checkpoint = torch.load(
    CHECKPOINT_PATH,
    map_location="cpu",
    weights_only=True
)

model.load_state_dict(
    checkpoint["model_state_dict"]
)

model.to(device)
model.eval()


# Last convolutional block.
target_layers = [
    model.layer4[-1]
]


transform = transforms.Compose([
    transforms.Resize(
        (224, 224)
    ),

    transforms.ToTensor(),

    transforms.Normalize(
        mean=[
            0.485,
            0.456,
            0.406
        ],

        std=[
            0.229,
            0.224,
            0.225
        ]
    )
])


# ============================================================
# Load paired analysis
# ============================================================

df = pd.read_csv(
    ERROR_PATH
)

df["id"] = (
    df["id"]
    .astype(str)
)


groups = [
    "fusion_only_correct",
    "roberta_only_correct",
    "both_correct",
    "both_wrong",
]


cam = GradCAM(
    model=model,
    target_layers=target_layers
)


summary_rows = []


for group in groups:

    subset = df[
        df["comparison_group"]
        == group
    ].copy()

    if len(subset) == 0:
        continue

    sample_n = min(
        N_PER_GROUP,
        len(subset)
    )

    sampled = subset.sample(
        n=sample_n,
        random_state=SEED
    )

    group_root = (
        OUTPUT_ROOT / group
    )

    group_root.mkdir(
        parents=True,
        exist_ok=True
    )


    print(
        "\n" + "=" * 70
    )

    print(
        group.upper()
    )

    print("=" * 70)


    for _, row in sampled.iterrows():

        image_path = Path(
            str(row["image_path"])
        )

        if not image_path.exists():

            print(
                "Missing:",
                image_path
            )

            continue


        with Image.open(
            image_path
        ) as image:

            image = image.convert(
                "RGB"
            )

            display_image = (
                image.resize(
                    (224, 224)
                )
            )

            rgb = (
                np.asarray(
                    display_image
                )
                .astype(np.float32)
                / 255.0
            )

            input_tensor = (
                transform(image)
                .unsqueeze(0)
                .to(device)
            )


        # Get ResNet's predicted class.
        with torch.no_grad():

            logits = model(
                input_tensor
            )

            predicted_class = int(
                torch.argmax(
                    logits,
                    dim=1
                ).item()
            )


        # Explain the predicted class.
        targets = [
            ClassifierOutputTarget(
                predicted_class
            )
        ]


        grayscale_cam = cam(
            input_tensor=input_tensor,
            targets=targets
        )[0]


        visualization = (
            show_cam_on_image(
                rgb,
                grayscale_cam,
                use_rgb=True
            )
        )


        output_path = (
            group_root
            / f"{row['id']}.jpg"
        )


        Image.fromarray(
            visualization
        ).save(
            output_path
        )


        summary_rows.append({
            "id":
                row["id"],

            "comparison_group":
                group,

            "label":
                int(row["label"]),

            "prediction_roberta":
                int(
                    row[
                        "prediction_roberta"
                    ]
                ),

            "prediction_resnet":
                int(
                    row[
                        "prediction_resnet"
                    ]
                ),

            "prediction_fusion":
                int(
                    row[
                        "prediction_fusion"
                    ]
                ),

            "probability_roberta":
                float(
                    row[
                        "probability_roberta"
                    ]
                ),

            "probability_resnet":
                float(
                    row[
                        "probability_resnet"
                    ]
                ),

            "probability_fused":
                float(
                    row[
                        "probability_fused"
                    ]
                ),

            "text":
                str(row["text"]),

            "image_path":
                str(image_path),

            "gradcam_path":
                str(output_path),
        })


        print(
            f"{row['id']} | "
            f"label={int(row['label'])} | "
            f"text={int(row['prediction_roberta'])} | "
            f"image={int(row['prediction_resnet'])} | "
            f"fusion={int(row['prediction_fusion'])}"
        )

# END REGISTERED SOURCE BLOCK


In [58]:
%%project_source multimodal-fake-news-detection/scripts/generate_gradcam_cases.py 1
summary = pd.DataFrame(
    summary_rows
)

summary.to_csv(
    OUTPUT_ROOT
    / "gradcam_case_summary.csv",
    index=False
)


print(
    "\n" + "=" * 70
)

print(
    "GRAD-CAM COMPLETE"
)

print("=" * 70)

print(
    f"\nGenerated {len(summary):,} "
    "case visualisations."
)

print(
    "Saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


### 6.7 Build multimodal case studies

Combine selected prediction and attribution evidence for inspection and reporting.

**Source:** `multimodal-fake-news-detection/scripts/build_multimodal_case_studies.py`  
**Imported modules:** `json`, `numpy`, `pandas`, `pathlib`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `results/gradcam/gradcam_case_summary.csv`
- `results/shap/all_token_attributions.csv`
- `results/case_studies`

The following cells contain the complete source; Run All registers it for inspection/export.

In [59]:
%%project_source multimodal-fake-news-detection/scripts/build_multimodal_case_studies.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd


GRADCAM_SUMMARY = Path(
    "results/gradcam/gradcam_case_summary.csv"
)

SHAP_TOKENS = Path(
    "results/shap/all_token_attributions.csv"
)

OUTPUT_ROOT = Path(
    "results/case_studies"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

N_PER_GROUP = 2

GROUPS = [
    "fusion_only_correct",
    "roberta_only_correct",
    "both_correct",
    "both_wrong",
]


# ============================================================
# Load Grad-CAM cases and SHAP token attributions
# ============================================================

gradcam = pd.read_csv(
    GRADCAM_SUMMARY
)

tokens = pd.read_csv(
    SHAP_TOKENS
)

gradcam["id"] = (
    gradcam["id"]
    .astype(str)
)

tokens["id"] = (
    tokens["id"]
    .astype(str)
)


# ============================================================
# Build corrected SHAP summaries
#
# Positive SHAP = supports explained RoBERTa class
# Negative SHAP = opposes explained RoBERTa class
# ============================================================

token_summaries = []


for sample_id, sample in tokens.groupby("id"):

        sample = sample[
        sample["token"].notna()
    ].copy()

        sample["token"] = (
        sample["token"]
        .astype(str)
    )

sample = sample[
        sample["token"]
        .str.strip()
        .ne("")
    ]


positive = (
        sample[
            sample["shap_value"] > 0
        ]
        .sort_values(
            "shap_value",
            ascending=False
        )
        .head(5)
    )

negative = (
        sample[
            sample["shap_value"] < 0
        ]
        .sort_values(
            "shap_value",
            ascending=True
        )
        .head(5)
    )


supportive = [
        {
            "token": str(row["token"]),
            "shap": float(
                row["shap_value"]
            ),
        }

        for _, row
        in positive.iterrows()
    ]


opposing = [
        {
            "token": str(row["token"]),
            "shap": float(
                row["shap_value"]
            ),
        }

        for _, row
        in negative.iterrows()
    ]


token_summaries.append({
        "id":
            sample_id,

        "supportive_tokens":
            json.dumps(
                supportive
            ),

        "opposing_tokens":
            json.dumps(
                opposing
            ),
    })


token_summary = pd.DataFrame(
    token_summaries
)


# ============================================================
# Merge SHAP + Grad-CAM case information
# ============================================================

df = gradcam.merge(
    token_summary,
    on="id",
    how="left",
    validate="one_to_one"
)


# ============================================================
# Calculate useful case-study characteristics
# ============================================================

# END REGISTERED SOURCE BLOCK


In [60]:
%%project_source multimodal-fake-news-detection/scripts/build_multimodal_case_studies.py 1
df["fusion_probability_shift"] = (
    df["probability_fused"]
    - df["probability_roberta"]
)

df["absolute_fusion_shift"] = (
    df["fusion_probability_shift"]
    .abs()
)


df["roberta_confidence"] = np.maximum(
    df["probability_roberta"],
    1.0 - df["probability_roberta"]
)

df["resnet_confidence"] = np.maximum(
    df["probability_resnet"],
    1.0 - df["probability_resnet"]
)

df["mean_model_confidence"] = (
    df["roberta_confidence"]
    + df["resnet_confidence"]
) / 2.0


# ============================================================
# Select two representative cases from each category
# ============================================================

selected_parts = []


for group in GROUPS:

    subset = df[
        df["comparison_group"]
        == group
    ].copy()


    if group in [
        "fusion_only_correct",
        "roberta_only_correct",
    ]:

        # For modality-conflict cases, select examples where
        # fusion moved the probability most strongly.
        subset = subset.sort_values(
            "absolute_fusion_shift",
            ascending=False
        )

    else:

        # For agreement / failure cases, select examples
        # where the unimodal models were most confident.
        subset = subset.sort_values(
            "mean_model_confidence",
            ascending=False
        )


    selected_parts.append(
        subset.head(
            N_PER_GROUP
        )
    )


selected = pd.concat(
    selected_parts,
    ignore_index=True
)


# ============================================================
# Save outputs
# ============================================================

df.to_csv(
    OUTPUT_ROOT
    / "all_32_multimodal_cases.csv",
    index=False
)

selected.to_csv(
    OUTPUT_ROOT
    / "selected_8_case_studies.csv",
    index=False
)


# ============================================================
# Print selected cases
# ============================================================

print("=" * 70)
print("MULTIMODAL CASE-STUDY CONSOLIDATION")
print("=" * 70)

print(
    f"\nAvailable explained cases: "
    f"{len(df)}"
)

print(
    f"Selected case studies: "
    f"{len(selected)}"
)


for group in GROUPS:

    group_df = selected[
        selected["comparison_group"]
        == group
    ]

    print(
        "\n" + "=" * 70
    )

    print(
        group.upper()
    )

    print("=" * 70)


    for _, row in group_df.iterrows():

        print(
            f"\nID: {row['id']}"
        )

        print(
            f"Text: {row['text']}"
        )

        print(
            f"True label: "
            f"{int(row['label'])}"
        )

        print(
            f"RoBERTa: "
            f"{int(row['prediction_roberta'])} "
            f"(P1={row['probability_roberta']:.3f})"
        )

        print(
            f"ResNet: "
            f"{int(row['prediction_resnet'])} "
            f"(P1={row['probability_resnet']:.3f})"
        )

        print(
            f"Fusion: "
            f"{int(row['prediction_fusion'])} "
            f"(P1={row['probability_fused']:.3f})"
        )

        print(
            "SHAP supporting:",
            row["supportive_tokens"]
        )

        print(
            "SHAP opposing:",
            row["opposing_tokens"]
        )

        print(
            "Grad-CAM:",
            row["gradcam_path"]
        )


# END REGISTERED SOURCE BLOCK


In [61]:
%%project_source multimodal-fake-news-detection/scripts/build_multimodal_case_studies.py 2
print(
    "\n" + "=" * 70
)

print(
    "CASE-STUDY CONSOLIDATION COMPLETE"
)

print("=" * 70)

print(
    "\nResults saved to:",
    OUTPUT_ROOT
)
# END REGISTERED SOURCE BLOCK


<a id="holdout"></a>
## 7. Locked final holdout

Do not repeatedly use this holdout to choose settings. Candidate construction, cleaning and freezing precede the final evaluation.

### 7.1 Create final holdout candidates

Select candidate cases for a separate final evaluation with the implemented exclusions.

**Source:** `multimodal-fake-news-detection/scripts/create_final_holdout_candidates.py`  
**Imported modules:** `json`, `pandas`, `pathlib`, `sklearn`  
**Top-level components:** `resolve_column`, `normalise_string`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/test.parquet`
- `data/processed/fakeddit/development`
- `data/processed/fakeddit/final_holdout`
- `results/metrics/final_holdout`

The following cells contain the complete source; Run All registers it for inspection/export.

In [62]:
%%project_source multimodal-fake-news-detection/scripts/create_final_holdout_candidates.py 0
import json
from pathlib import Path

import pandas as pd
from sklearn.model_selection import train_test_split


SEED = 2026
CANDIDATE_SIZE = 10000


FULL_TEST_PATH = Path(
    "data/processed/fakeddit/test.parquet"
)

DEV_ROOT = Path(
    "data/processed/fakeddit/development"
)

OUTPUT_ROOT = Path(
    "data/processed/fakeddit/final_holdout"
)

METRICS_ROOT = Path(
    "results/metrics/final_holdout"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

METRICS_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


def resolve_column(
    dataframe,
    candidates,
    name
):

    for column in candidates:

        if column in dataframe.columns:
            return column

    raise ValueError(
        f"Could not find {name}. "
        f"Available columns: "
        f"{list(dataframe.columns)}"
    )


def normalise_string(series):

    return (
        series
        .astype("string")
        .fillna("")
        .str.strip()
    )


print("=" * 70)
print("CREATE FINAL HOLDOUT CANDIDATES")
print("=" * 70)


# ============================================================
# Load full official public test pool
# ============================================================

full = pd.read_parquet(
    FULL_TEST_PATH
)

print(
    f"\nFull public test rows: "
    f"{len(full):,}"
)

print(
    "\nColumns:"
)

print(
    list(full.columns)
)


id_col = resolve_column(
    full,
    ["id"],
    "ID column"
)

label_col = resolve_column(
    full,
    [
        "label",
        "2_way_label",
    ],
    "binary label column"
)

text_col = resolve_column(
    full,
    [
        "text",
        "clean_title",
        "title",
    ],
    "text column"
)

image_url_col = resolve_column(
    full,
    [
        "image_url",
    ],
    "image URL column"
)


# ============================================================
# Load ALL development manifests
#
# These include every sample we have previously used:
# train + validation + development test.
# ============================================================

development_frames = []

for split in [
    "train",
    "validation",
    "test",
]:

    path = (
        DEV_ROOT
        / f"{split}.parquet"
    )

    frame = pd.read_parquet(
        path
    )

    frame["_development_split"] = (
        split
    )

    development_frames.append(
        frame
    )


# END REGISTERED SOURCE BLOCK


In [63]:
%%project_source multimodal-fake-news-detection/scripts/create_final_holdout_candidates.py 1
development = pd.concat(
    development_frames,
    ignore_index=True
)


print(
    f"\nPreviously used development rows: "
    f"{len(development):,}"
)


dev_id_col = resolve_column(
    development,
    ["id"],
    "development ID column"
)

dev_text_col = resolve_column(
    development,
    [
        "text",
        "clean_title",
        "title",
    ],
    "development text column"
)

dev_image_url_col = resolve_column(
    development,
    ["image_url"],
    "development image URL column"
)


# ============================================================
# Canonical values for overlap checks
# ============================================================

full_ids = normalise_string(
    full[id_col]
)

full_text = normalise_string(
    full[text_col]
)

full_urls = normalise_string(
    full[image_url_col]
)


development_ids = set(
    normalise_string(
        development[dev_id_col]
    )
)

development_text = set(
    value
    for value in normalise_string(
        development[dev_text_col]
    )
    if value != ""
)

development_urls = set(
    value
    for value in normalise_string(
        development[dev_image_url_col]
    )
    if value != ""
)


# ============================================================
# Leakage exclusion
#
# Final holdout cannot share:
# - ID
# - exact processed text
# - exact image URL
#
# with anything previously used during development.
# ============================================================

id_overlap = (
    full_ids.isin(
        development_ids
    )
)

text_overlap = (
    full_text.ne("")
    &
    full_text.isin(
        development_text
    )
)

url_overlap = (
    full_urls.ne("")
    &
    full_urls.isin(
        development_urls
    )
)


any_overlap = (
    id_overlap
    |
    text_overlap
    |
    url_overlap
)


print(
    "\nOverlap with development data:"
)

print(
    f"ID overlap:        "
    f"{int(id_overlap.sum()):,}"
)

print(
    f"Exact text overlap:"
    f" {int(text_overlap.sum()):,}"
)

print(
    f"Image URL overlap: "
    f"{int(url_overlap.sum()):,}"
)

print(
    f"Excluded by union: "
    f"{int(any_overlap.sum()):,}"
)


eligible = (
    full.loc[
        ~any_overlap
    ]
    .copy()
    .reset_index(drop=True)
)


print(
    f"\nEligible untouched pool: "
    f"{len(eligible):,}"
)


if len(eligible) < CANDIDATE_SIZE:

    raise ValueError(
        "Eligible pool is smaller than "
        f"{CANDIDATE_SIZE:,}."
    )


# ============================================================
# Select 10,000 candidates
#
# Stratification preserves the binary-label distribution
# of the untouched eligible pool.
# ============================================================

# END REGISTERED SOURCE BLOCK


In [64]:
%%project_source multimodal-fake-news-detection/scripts/create_final_holdout_candidates.py 2
candidates, _ = train_test_split(
    eligible,
    train_size=CANDIDATE_SIZE,
    random_state=SEED,
    stratify=eligible[label_col],
)


candidates = (
    candidates
    .sample(
        frac=1.0,
        random_state=SEED
    )
    .reset_index(drop=True)
)


# Standard aliases for downstream scripts.
candidates["id"] = (
    candidates[id_col]
    .astype(str)
)

candidates["label"] = (
    candidates[label_col]
    .astype(int)
)

candidates["text"] = (
    candidates[text_col]
    .astype("string")
    .fillna("")
)

candidates["image_url"] = (
    candidates[image_url_col]
    .astype("string")
    .fillna("")
)


output_path = (
    OUTPUT_ROOT
    / "candidates.parquet"
)

candidates.to_parquet(
    output_path,
    index=False
)


# ============================================================
# Reproducibility metadata
# ============================================================

label_counts = {
    str(key): int(value)
    for key, value
    in candidates[
        "label"
    ]
    .value_counts()
    .sort_index()
    .items()
}


metadata = {
    "purpose":
        "unseen final evaluation holdout",

    "source":
        str(FULL_TEST_PATH),

    "candidate_seed":
        SEED,

    "candidate_size":
        CANDIDATE_SIZE,

    "full_public_test_rows":
        int(len(full)),

    "previous_development_rows":
        int(len(development)),

    "overlap_counts": {
        "id":
            int(id_overlap.sum()),

        "exact_text":
            int(text_overlap.sum()),

        "image_url":
            int(url_overlap.sum()),

        "union_excluded":
            int(any_overlap.sum()),
    },

    "eligible_pool_rows":
        int(len(eligible)),

    "candidate_label_counts":
        label_counts,

    "model_predictions_used":
        False,

    "test_metrics_used_for_selection":
        False,
}


with (
    METRICS_ROOT
    / "candidate_selection.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        metadata,
        f,
        indent=2
    )


print(
    "\nCandidate label counts:"
)

print(
    candidates[
        "label"
    ]
    .value_counts()
    .sort_index()
)


print(
    "\nCandidate manifest saved to:"
)

print(
    output_path
)


print(
    "\nIMPORTANT:"
)

print(
    "No model predictions or model "
    "performance were used to select "
    "these samples."
)


# END REGISTERED SOURCE BLOCK


In [65]:
%%project_source multimodal-fake-news-detection/scripts/create_final_holdout_candidates.py 3
print(
    "\n" + "=" * 70
)

print(
    "FINAL HOLDOUT CANDIDATE "
    "SELECTION COMPLETE"
)

print("=" * 70)
# END REGISTERED SOURCE BLOCK


### 7.2 Prepare final holdout

Acquire and audit final candidate images, exclude invalid content and prepare the locked usable holdout records.

**Source:** `multimodal-fake-news-detection/scripts/prepare_final_holdout.py`  
**Imported modules:** `PIL`, `concurrent`, `hashlib`, `io`, `json`, `pandas`, `pathlib`, `requests`, `time`  
**Top-level components:** `sha256_bytes`, `sha256_file`, `validate_image_bytes`, `validate_existing_file`, `download_one`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/final_holdout/candidates.parquet`
- `data/raw/fakeddit/final_holdout_images`
- `data/raw/fakeddit/development_images`
- `data/processed/fakeddit/final_holdout`
- `results/metrics/final_holdout`

The following cells contain the complete source; Run All registers it for inspection/export.

In [66]:
%%project_source multimodal-fake-news-detection/scripts/prepare_final_holdout.py 0
import hashlib
import json
import time
from concurrent.futures import ThreadPoolExecutor, as_completed
from io import BytesIO
from pathlib import Path

import pandas as pd
import requests
from PIL import Image


CANDIDATE_PATH = Path(
    "data/processed/fakeddit/final_holdout/candidates.parquet"
)

IMAGE_ROOT = Path(
    "data/raw/fakeddit/final_holdout_images"
)

DEVELOPMENT_IMAGE_ROOT = Path(
    "data/raw/fakeddit/development_images"
)

OUTPUT_ROOT = Path(
    "data/processed/fakeddit/final_holdout"
)

METRICS_ROOT = Path(
    "results/metrics/final_holdout"
)


FINAL_SIZE = 5000

MAX_WORKERS = 16
TIMEOUT_SECONDS = 20
MAX_ATTEMPTS = 3


# Known invalid "not available in your region" placeholder.
PLACEHOLDER_HASH = (
    "faa24ec881e6040655c187a681d6dc496eb8aa41e1bd0652a180b3a40b457187"
)


IMAGE_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)

METRICS_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


HEADERS = {
    "User-Agent":
        "Mozilla/5.0 multimodal-fake-news-research"
}


def sha256_bytes(data):

    return hashlib.sha256(
        data
    ).hexdigest()


def sha256_file(path):

    digest = hashlib.sha256()

    with path.open("rb") as f:

        for chunk in iter(
            lambda: f.read(1024 * 1024),
            b""
        ):
            digest.update(chunk)

    return digest.hexdigest()


def validate_image_bytes(data):

    try:

        with Image.open(
            BytesIO(data)
        ) as image:

            image.verify()

        # Open a second time because verify()
        # invalidates the first PIL object.
        with Image.open(
            BytesIO(data)
        ) as image:

            image = image.convert("RGB")

            width, height = image.size

        return (
            True,
            int(width),
            int(height),
            None,
        )

    except Exception as exc:

        return (
            False,
            None,
            None,
            str(exc),
        )


def validate_existing_file(path):

    try:

        data = path.read_bytes()

    except Exception as exc:

        return {
            "valid":
                False,

            "sha256":
                None,

            "width":
                None,

            "height":
                None,

            "error":
                str(exc),
        }


    valid, width, height, error = (
        validate_image_bytes(data)
    )

    return {
        "valid":
            valid,

        "sha256":
            (
                sha256_bytes(data)
                if valid
                else None
            ),

        "width":
            width,

        "height":
            height,

        "error":
            error,
    }


# END REGISTERED SOURCE BLOCK


In [67]:
%%project_source multimodal-fake-news-detection/scripts/prepare_final_holdout.py 1
def download_one(index, row):

    sample_id = str(
        row["id"]
    )

    url = str(
        row["image_url"]
    ).strip()

    output_path = (
        IMAGE_ROOT
        / f"{sample_id}.jpg"
    )


    result = {
        "candidate_order":
            int(index),

        "id":
            sample_id,

        "image_path":
            str(output_path),

        "download_status":
            None,

        "image_valid":
            False,

        "image_sha256":
            None,

        "image_width":
            None,

        "image_height":
            None,

        "download_error":
            None,
    }


    if (
        not url
        or url.lower() == "nan"
    ):

        result[
            "download_status"
        ] = "missing_url"

        return result


    # --------------------------------------------------------
    # Reuse an existing downloaded file.
    # --------------------------------------------------------

    if output_path.exists():

        checked = (
            validate_existing_file(
                output_path
            )
        )

        if checked["valid"]:

            result.update({
                "download_status":
                    "already_present",

                "image_valid":
                    True,

                "image_sha256":
                    checked["sha256"],

                "image_width":
                    checked["width"],

                "image_height":
                    checked["height"],
            })

            return result

        else:

            # Remove broken partial download
            # and try again.
            try:
                output_path.unlink()
            except Exception:
                pass


    # --------------------------------------------------------
    # Download with retry.
    # --------------------------------------------------------

    last_error = None


    for attempt in range(
        1,
        MAX_ATTEMPTS + 1
    ):

        try:

            response = requests.get(
                url,
                headers=HEADERS,
                timeout=TIMEOUT_SECONDS
            )

            response.raise_for_status()

            data = response.content


            valid, width, height, error = (
                validate_image_bytes(
                    data
                )
            )


            if not valid:

                last_error = (
                    f"invalid_image: {error}"
                )

                continue


            output_path.write_bytes(
                data
            )


            result.update({
                "download_status":
                    "downloaded",

                "image_valid":
                    True,

                "image_sha256":
                    sha256_bytes(data),

                "image_width":
                    width,

                "image_height":
                    height,

                "download_error":
                    None,
            })


            return result


        except Exception as exc:

            last_error = str(exc)

            if attempt < MAX_ATTEMPTS:

                time.sleep(
                    0.5 * attempt
                )


    result[
        "download_status"
    ] = "failed"

    result[
        "download_error"
    ] = last_error

    return result


# END REGISTERED SOURCE BLOCK


In [68]:
%%project_source multimodal-fake-news-detection/scripts/prepare_final_holdout.py 2
print("=" * 70)
print("PREPARE FINAL UNSEEN HOLDOUT")
print("=" * 70)


# ============================================================
# Load frozen candidate manifest
# ============================================================

candidates = pd.read_parquet(
    CANDIDATE_PATH
)

candidates["id"] = (
    candidates["id"]
    .astype(str)
)

candidates["text"] = (
    candidates["text"]
    .astype("string")
    .fillna("")
)

candidates["image_url"] = (
    candidates["image_url"]
    .astype("string")
    .fillna("")
)


print(
    f"\nFrozen candidates: "
    f"{len(candidates):,}"
)

print(
    f"Target final holdout: "
    f"{FINAL_SIZE:,}"
)


# ============================================================
# Hash all EXISTING development images
#
# This detects visual duplicates even when URLs differ.
# ============================================================

print(
    "\nHashing existing development images..."
)


development_hashes = set()

development_files = [
    path
    for path
    in DEVELOPMENT_IMAGE_ROOT.rglob("*")
    if path.is_file()
]


for i, path in enumerate(
    development_files,
    start=1
):

    try:

        development_hashes.add(
            sha256_file(path)
        )

    except Exception:
        pass


    if i % 5000 == 0:

        print(
            f"  Hashed {i:,} "
            "development files"
        )


print(
    f"Development files scanned: "
    f"{len(development_files):,}"
)

print(
    f"Unique development image hashes: "
    f"{len(development_hashes):,}"
)


# ============================================================
# Download candidate images
# ============================================================

print(
    "\nDownloading / validating "
    "candidate images..."
)

print(
    f"Workers: {MAX_WORKERS}"
)


records = []


with ThreadPoolExecutor(
    max_workers=MAX_WORKERS
) as executor:

    futures = {
        executor.submit(
            download_one,
            index,
            row
        ): index

        for index, row
        in candidates.iterrows()
    }


    completed = 0


    for future in as_completed(
        futures
    ):

        records.append(
            future.result()
        )

        completed += 1


        if (
            completed % 500 == 0
            or completed
            == len(candidates)
        ):

            print(
                f"  Completed "
                f"{completed:,} / "
                f"{len(candidates):,}"
            )


status = pd.DataFrame(
    records
)


# Restore deterministic candidate order.
# END REGISTERED SOURCE BLOCK


In [69]:
%%project_source multimodal-fake-news-detection/scripts/prepare_final_holdout.py 3
status = status.sort_values(
    "candidate_order"
).reset_index(
    drop=True
)


manifest = candidates.merge(
    status,
    on="id",
    how="left",
    validate="one_to_one"
)


# ============================================================
# Cleaning flags
# ============================================================

manifest[
    "is_known_placeholder"
] = (
    manifest["image_sha256"]
    == PLACEHOLDER_HASH
)


manifest[
    "image_seen_in_development"
] = (
    manifest["image_sha256"]
    .fillna("")
    .isin(
        development_hashes
    )
)


# Exact duplicate text within final candidate pool.
#
# Keep the earliest sample in the already-frozen
# candidate order.
normalised_text = (
    manifest["text"]
    .astype("string")
    .fillna("")
    .str.strip()
)

manifest[
    "duplicate_text_within_candidates"
] = (
    normalised_text.ne("")
    &
    normalised_text.duplicated(
        keep="first"
    )
)


# Exact image duplicate inside final candidate pool.
#
# Again keep first occurrence only.
hash_values = (
    manifest[
        "image_sha256"
    ]
    .fillna("")
)

manifest[
    "duplicate_image_within_candidates"
] = (
    hash_values.ne("")
    &
    hash_values.duplicated(
        keep="first"
    )
)


manifest[
    "usable_final"
] = (
    manifest[
        "image_valid"
    ].fillna(False)
    &
    ~manifest[
        "is_known_placeholder"
    ]
    &
    ~manifest[
        "image_seen_in_development"
    ]
    &
    ~manifest[
        "duplicate_text_within_candidates"
    ]
    &
    ~manifest[
        "duplicate_image_within_candidates"
    ]
)


# ============================================================
# Diagnostics
# ============================================================

print(
    "\nDownload status:"
)

print(
    manifest[
        "download_status"
    ]
    .value_counts(
        dropna=False
    )
)


print(
    "\nCleaning exclusions:"
)

print(
    "Invalid / unavailable image:",
    int(
        (
            ~manifest[
                "image_valid"
            ].fillna(False)
        ).sum()
    )
)

print(
    "Known placeholder:",
    int(
        manifest[
            "is_known_placeholder"
        ].sum()
    )
)

print(
    "Image seen in development:",
    int(
        manifest[
            "image_seen_in_development"
        ].sum()
    )
)

print(
    "Duplicate text within candidates:",
    int(
        manifest[
            "duplicate_text_within_candidates"
        ].sum()
    )
)

# END REGISTERED SOURCE BLOCK


In [70]:
%%project_source multimodal-fake-news-detection/scripts/prepare_final_holdout.py 4
print(
    "Duplicate image within candidates:",
    int(
        manifest[
            "duplicate_image_within_candidates"
        ].sum()
    )
)


usable = manifest[
    manifest[
        "usable_final"
    ]
].copy()


print(
    f"\nUsable leakage-reduced samples: "
    f"{len(usable):,}"
)


if len(usable) < FINAL_SIZE:

    raise RuntimeError(
        "Fewer than "
        f"{FINAL_SIZE:,} usable samples. "
        "Do not change model settings. "
        "Increase the candidate pool instead."
    )


# ============================================================
# Freeze EXACTLY first 5,000 usable samples
#
# Candidate ordering was fixed before any image download
# or model evaluation.
# ============================================================

final = (
    usable
    .head(
        FINAL_SIZE
    )
    .copy()
    .reset_index(drop=True)
)


# ============================================================
# Final overlap assertions
# ============================================================

assert (
    final["id"]
    .nunique()
    == len(final)
)

assert not final[
    "is_known_placeholder"
].any()

assert not final[
    "image_seen_in_development"
].any()

assert not final[
    "duplicate_text_within_candidates"
].any()

assert not final[
    "duplicate_image_within_candidates"
].any()


# ============================================================
# Holdout fingerprint
# ============================================================

ordered_ids = "\n".join(
    final["id"]
    .astype(str)
    .tolist()
)

id_sha256 = hashlib.sha256(
    ordered_ids.encode("utf-8")
).hexdigest()


# ============================================================
# Save manifests
# ============================================================

manifest.to_parquet(
    OUTPUT_ROOT
    / "candidate_image_status.parquet",
    index=False
)

final.to_parquet(
    OUTPUT_ROOT
    / "final_5000.parquet",
    index=False
)


label_counts = {
    str(key): int(value)
    for key, value
    in final[
        "label"
    ]
    .value_counts()
    .sort_index()
    .items()
}


metadata = {
    "purpose":
        "final unseen multimodal evaluation",

    "candidate_count":
        int(len(candidates)),

    "target_final_count":
        FINAL_SIZE,

    "usable_before_final_selection":
        int(len(usable)),

    "final_count":
        int(len(final)),

    "final_label_counts":
        label_counts,

    "ordered_id_sha256":
        id_sha256,

    "known_placeholder_hash":
        PLACEHOLDER_HASH,

    "cleaning": {
        "require_readable_image":
            True,

        "exclude_known_placeholder":
            True,

        "exclude_development_image_hashes":
            True,

        "deduplicate_exact_text_within_candidates":
            True,

        "deduplicate_exact_image_hash_within_candidates":
            True,
    },

    "fusion_model_locked": {
        "text_model":
            "roberta-base fine-tuned checkpoint",

        "image_model":
            "resnet50 fine-tuned checkpoint",

        "alpha_text":
            0.45,

        "alpha_image":
            0.55,

        "decision_threshold":
            0.5,
    },

    "model_predictions_used_for_selection":
        False,

    "model_metrics_used_for_selection":
        False,
}


# END REGISTERED SOURCE BLOCK


In [71]:
%%project_source multimodal-fake-news-detection/scripts/prepare_final_holdout.py 5
with (
    METRICS_ROOT
    / "final_holdout_freeze.json"
).open(
    "w",
    encoding="utf-8"
) as f:

    json.dump(
        metadata,
        f,
        indent=2
    )


print(
    "\n" + "=" * 70
)

print(
    "FINAL HOLDOUT FROZEN"
)

print("=" * 70)


print(
    f"\nFinal samples: "
    f"{len(final):,}"
)

print(
    "\nFinal label counts:"
)

print(
    final[
        "label"
    ]
    .value_counts()
    .sort_index()
)


print(
    "\nOrdered ID SHA256:"
)

print(
    id_sha256
)


print(
    "\nFinal manifest:"
)

print(
    OUTPUT_ROOT
    / "final_5000.parquet"
)


print(
    "\nIMPORTANT:"
)

print(
    "The final holdout is now frozen."
)

print(
    "Do not alter models, fusion weights, "
    "thresholds, or cleaning rules after "
    "viewing final performance."
)
# END REGISTERED SOURCE BLOCK


### 7.3 Evaluate final holdout

Apply frozen settings to the final holdout, record predictions, metrics, paired comparisons and calibration.

**Source:** `multimodal-fake-news-detection/scripts/evaluate_final_holdout.py`  
**Imported modules:** `PIL`, `hashlib`, `json`, `numpy`, `pandas`, `pathlib`, `scipy`, `sklearn`, `torch`, `torchvision`, `transformers`  
**Top-level components:** `TextDataset`, `ImageDataset`, `calculate_metrics`, `expected_calibration_error`, `predict_roberta`, `predict_resnet`, `paired_bootstrap`, `main`

**Literal data/output path references** (inspect the code for read/write direction and constructed paths):
- `data/processed/fakeddit/final_holdout/final_5000.parquet`
- `checkpoints/roberta_baseline`
- `checkpoints/resnet50_baseline/best_model.pt`
- `results/metrics/final_evaluation`

The following cells contain the complete source; Run All registers it for inspection/export.

In [72]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_final_holdout.py 0
import json
from pathlib import Path

import numpy as np
import pandas as pd
from PIL import Image

import torch
import torch.nn as nn
from torch.utils.data import Dataset, DataLoader

from transformers import (
    AutoTokenizer,
    AutoModelForSequenceClassification,
)

from torchvision.models import resnet50
from torchvision import transforms

from sklearn.metrics import (
    accuracy_score,
    precision_score,
    recall_score,
    f1_score,
    roc_auc_score,
    average_precision_score,
    confusion_matrix,
    brier_score_loss,
    log_loss,
)

from scipy.stats import binomtest


# ============================================================
# LOCKED FINAL SPECIFICATION
# ============================================================

FINAL_MANIFEST = Path(
    "data/processed/fakeddit/final_holdout/final_5000.parquet"
)

ROBERTA_CHECKPOINT = Path(
    "checkpoints/roberta_baseline"
)

RESNET_CHECKPOINT = Path(
    "checkpoints/resnet50_baseline/best_model.pt"
)

OUTPUT_ROOT = Path(
    "results/metrics/final_evaluation"
)

OUTPUT_ROOT.mkdir(
    parents=True,
    exist_ok=True
)


ALPHA_TEXT = 0.45
ALPHA_IMAGE = 0.55

THRESHOLD = 0.50

MAX_LENGTH = 64

ROBERTA_BATCH_SIZE = 16
RESNET_BATCH_SIZE = 32

NUM_WORKERS = 4

BOOTSTRAP_SAMPLES = 5000
BOOTSTRAP_SEED = 42

EXPECTED_HOLDOUT_SIZE = 5000

EXPECTED_ID_SHA256 = (
    "2ebe8ee8bf208f291f65c67c069e38a2922ec89af80387d94a865417a914494a"
)


# ============================================================
# Dataset classes
# ============================================================

class TextDataset(Dataset):

    def __init__(
        self,
        dataframe,
        tokenizer
    ):

        self.df = (
            dataframe
            .reset_index(drop=True)
        )

        self.tokenizer = tokenizer


    def __len__(self):

        return len(self.df)


    def __getitem__(
        self,
        idx
    ):

        row = self.df.iloc[idx]

        encoded = self.tokenizer(
            str(row["text"]),
            padding="max_length",
            truncation=True,
            max_length=MAX_LENGTH,
            return_tensors="pt"
        )

        return {
            "id":
                str(row["id"]),

            "label":
                int(row["label"]),

            "input_ids":
                encoded[
                    "input_ids"
                ].squeeze(0),

            "attention_mask":
                encoded[
                    "attention_mask"
                ].squeeze(0),
        }


class ImageDataset(Dataset):

    def __init__(
        self,
        dataframe,
        transform
    ):

        self.df = (
            dataframe
            .reset_index(drop=True)
        )

        self.transform = transform


    def __len__(self):

        return len(self.df)


    def __getitem__(
        self,
        idx
    ):

        row = self.df.iloc[idx]

        image_path = Path(
            str(row["image_path"])
        )

        with Image.open(
            image_path
        ) as image:

            image = image.convert(
                "RGB"
            )

            image = self.transform(
                image
            )

        return {
            "id":
                str(row["id"]),

            "label":
                int(row["label"]),

            "image":
                image,
        }


# ============================================================
# Metrics
# ============================================================

# END REGISTERED SOURCE BLOCK


In [73]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_final_holdout.py 1
def calculate_metrics(
    labels,
    predictions,
    probabilities
):

    return {
        "accuracy":
            float(
                accuracy_score(
                    labels,
                    predictions
                )
            ),

        "precision":
            float(
                precision_score(
                    labels,
                    predictions,
                    zero_division=0
                )
            ),

        "recall":
            float(
                recall_score(
                    labels,
                    predictions,
                    zero_division=0
                )
            ),

        "f1":
            float(
                f1_score(
                    labels,
                    predictions,
                    zero_division=0
                )
            ),

        "f1_macro":
            float(
                f1_score(
                    labels,
                    predictions,
                    average="macro",
                    zero_division=0
                )
            ),

        "roc_auc":
            float(
                roc_auc_score(
                    labels,
                    probabilities
                )
            ),

        "pr_auc":
            float(
                average_precision_score(
                    labels,
                    probabilities
                )
            ),

        "brier_score":
            float(
                brier_score_loss(
                    labels,
                    probabilities
                )
            ),

        "log_loss":
            float(
                log_loss(
                    labels,
                    np.clip(
                        probabilities,
                        1e-7,
                        1 - 1e-7
                    )
                )
            ),

        "confusion_matrix":
            confusion_matrix(
                labels,
                predictions
            ).tolist(),
    }


def expected_calibration_error(
    labels,
    probabilities,
    n_bins=10
):

    labels = np.asarray(
        labels
    )

    probabilities = np.asarray(
        probabilities
    )

    predictions = (
        probabilities
        >= THRESHOLD
    ).astype(int)

    confidence = np.maximum(
        probabilities,
        1.0 - probabilities
    )

    correctness = (
        predictions
        == labels
    ).astype(float)

    edges = np.linspace(
        0.5,
        1.0,
        n_bins + 1
    )

    ece = 0.0


    for i in range(
        n_bins
    ):

        lower = edges[i]
        upper = edges[i + 1]

        if i == n_bins - 1:

            mask = (
                (confidence >= lower)
                &
                (confidence <= upper)
            )

        else:

            mask = (
                (confidence >= lower)
                &
                (confidence < upper)
            )


        if not mask.any():
            continue


        bin_accuracy = (
            correctness[
                mask
            ].mean()
        )

        bin_confidence = (
            confidence[
                mask
            ].mean()
        )


        ece += (
            mask.mean()
            *
            abs(
                bin_accuracy
                - bin_confidence
            )
        )


    return float(ece)


# ============================================================
# Inference
# ============================================================

# END REGISTERED SOURCE BLOCK


In [74]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_final_holdout.py 2
@torch.no_grad()
def predict_roberta(
    dataframe,
    model,
    tokenizer,
    device
):

    dataset = TextDataset(
        dataframe,
        tokenizer
    )

    loader = DataLoader(
        dataset,
        batch_size=ROBERTA_BATCH_SIZE,
        shuffle=False,
        num_workers=0,
        pin_memory=(
            device.type
            == "cuda"
        )
    )

    ids = []
    labels = []
    probabilities = []


    model.eval()


    for batch in loader:

        input_ids = (
            batch[
                "input_ids"
            ]
            .to(
                device,
                non_blocking=True
            )
        )

        attention_mask = (
            batch[
                "attention_mask"
            ]
            .to(
                device,
                non_blocking=True
            )
        )


        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=(
                device.type
                == "cuda"
            )
        ):

            logits = model(
                input_ids=input_ids,
                attention_mask=attention_mask
            ).logits


        probs = torch.softmax(
            logits,
            dim=1
        )[:, 1]


        ids.extend(
            batch["id"]
        )

        labels.extend(
            batch["label"]
            .numpy()
            .tolist()
        )

        probabilities.extend(
            probs
            .cpu()
            .numpy()
            .tolist()
        )


    probabilities = np.asarray(
        probabilities
    )

    predictions = (
        probabilities
        >= THRESHOLD
    ).astype(int)


    return pd.DataFrame({
        "id":
            ids,

        "label":
            labels,

        "probability_roberta":
            probabilities,

        "prediction_roberta":
            predictions,
    })


@torch.no_grad()
def predict_resnet(
    dataframe,
    model,
    transform,
    device
):

    dataset = ImageDataset(
        dataframe,
        transform
    )


    loader_kwargs = {
        "batch_size":
            RESNET_BATCH_SIZE,

        "shuffle":
            False,

        "num_workers":
            NUM_WORKERS,

        "pin_memory":
            (
                device.type
                == "cuda"
            ),
    }


    if NUM_WORKERS > 0:

        loader_kwargs[
            "persistent_workers"
        ] = True


    loader = DataLoader(
        dataset,
        **loader_kwargs
    )


    ids = []
    labels = []
    probabilities = []


    model.eval()


    for batch in loader:

        images = (
            batch["image"]
            .to(
                device,
                non_blocking=True
            )
        )


        with torch.autocast(
            device_type="cuda",
            dtype=torch.float16,
            enabled=(
                device.type
                == "cuda"
            )
        ):

            logits = model(
                images
            )


        probs = torch.softmax(
            logits,
            dim=1
        )[:, 1]


        ids.extend(
            batch["id"]
        )

        labels.extend(
            batch["label"]
            .numpy()
            .tolist()
        )

        probabilities.extend(
            probs
            .cpu()
            .numpy()
            .tolist()
        )


    probabilities = np.asarray(
        probabilities
    )

    predictions = (
        probabilities
        >= THRESHOLD
    ).astype(int)


    return pd.DataFrame({
        "id":
            ids,

        "label":
            labels,

        "probability_resnet":
            probabilities,

        "prediction_resnet":
            predictions,
    })


# ============================================================
# Paired bootstrap
# ============================================================

# END REGISTERED SOURCE BLOCK


In [75]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_final_holdout.py 3
def paired_bootstrap(
    labels,
    baseline_pred,
    baseline_prob,
    fusion_pred,
    fusion_prob
):

    rng = np.random.default_rng(
        BOOTSTRAP_SEED
    )

    n = len(labels)


    metric_names = [
        "accuracy",
        "f1",
        "f1_macro",
        "roc_auc",
        "pr_auc",
    ]


    differences = {
        metric: []
        for metric
        in metric_names
    }


    for _ in range(
        BOOTSTRAP_SAMPLES
    ):

        indices = rng.integers(
            0,
            n,
            size=n
        )

        y_sample = labels[
            indices
        ]


        if (
            len(
                np.unique(
                    y_sample
                )
            )
            < 2
        ):
            continue


        baseline = calculate_metrics(
            y_sample,
            baseline_pred[
                indices
            ],
            baseline_prob[
                indices
            ]
        )

        fused = calculate_metrics(
            y_sample,
            fusion_pred[
                indices
            ],
            fusion_prob[
                indices
            ]
        )


        for metric in metric_names:

            differences[
                metric
            ].append(
                fused[metric]
                -
                baseline[metric]
            )


    output = {}


    for metric in metric_names:

        values = np.asarray(
            differences[
                metric
            ]
        )

        output[
            metric
        ] = {
            "ci_95_lower":
                float(
                    np.percentile(
                        values,
                        2.5
                    )
                ),

            "ci_95_upper":
                float(
                    np.percentile(
                        values,
                        97.5
                    )
                ),
        }


    return output


# ============================================================
# Main
# ============================================================

def main():

    print("=" * 70)
    print("FINAL UNSEEN HOLDOUT EVALUATION")
    print("=" * 70)


    dataframe = pd.read_parquet(
        FINAL_MANIFEST
    )


    if (
        len(dataframe)
        != EXPECTED_HOLDOUT_SIZE
    ):

        raise ValueError(
            "Final holdout size mismatch."
        )


    # Verify exact ordered holdout fingerprint.
    import hashlib

    ordered_ids = "\n".join(
        dataframe[
            "id"
        ]
        .astype(str)
        .tolist()
    )

    fingerprint = hashlib.sha256(
        ordered_ids.encode(
            "utf-8"
        )
    ).hexdigest()


    print(
        f"\nSamples: "
        f"{len(dataframe):,}"
    )

    print(
        "Holdout SHA256:",
        fingerprint
    )


    if (
        fingerprint
        != EXPECTED_ID_SHA256
    ):

        raise ValueError(
            "FINAL HOLDOUT FINGERPRINT "
            "DOES NOT MATCH LOCKED SET."
        )


    print(
        "\nHoldout fingerprint verified."
    )


    print(
        "\nLabel counts:"
    )

    print(
        dataframe[
            "label"
        ]
        .value_counts()
        .sort_index()
    )


    device = torch.device(
        "cuda"
        if torch.cuda.is_available()
        else "cpu"
    )


    print(
        f"\nDevice: {device}"
    )

    if (
        device.type
        == "cuda"
    ):

        print(
            "GPU:",
            torch.cuda.get_device_name(
                0
            )
        )


    # ========================================================
    # Load locked RoBERTa
    # ========================================================

    print(
        "\nLoading locked RoBERTa..."
    )

    tokenizer = (
        AutoTokenizer
        .from_pretrained(
            ROBERTA_CHECKPOINT
        )
    )

    roberta = (
        AutoModelForSequenceClassification
        .from_pretrained(
            ROBERTA_CHECKPOINT
        )
    )

    roberta.to(
        device
    )


    # ========================================================
    # Load locked ResNet
    # ========================================================

    print(
        "Loading locked ResNet..."
    )

    checkpoint = torch.load(
        RESNET_CHECKPOINT,
        map_location="cpu",
        weights_only=True
    )

    resnet = resnet50(
        weights=None
    )

    features = (
        resnet.fc.in_features
    )

    resnet.fc = nn.Linear(
        features,
        2
    )

    resnet.load_state_dict(
        checkpoint[
            "model_state_dict"
        ]
    )

    resnet.to(
        device
    )


    image_transform = transforms.Compose([
        transforms.Resize(
            (224, 224)
        ),

        transforms.ToTensor(),

        transforms.Normalize(
            mean=[
                0.485,
                0.456,
                0.406,
            ],

            std=[
                0.229,
                0.224,
                0.225,
            ]
        ),
    ])


    # ========================================================
    # FINAL inference
    # ========================================================

    print(
        "\nRunning RoBERTa inference..."
    )

    text_results = predict_roberta(
        dataframe,
        roberta,
        tokenizer,
        device
    )


    print(
        "Running ResNet inference..."
    )

    image_results = predict_resnet(
        dataframe,
        resnet,
        image_transform,
        device
    )


    results = text_results.merge(
        image_results[
            [
                "id",
                "probability_resnet",
                "prediction_resnet",
            ]
        ],
        on="id",
        validate="one_to_one"
    )


    # ========================================================
    # LOCKED late fusion
    # ========================================================

    results[
        "probability_fusion"
    ] = (
        ALPHA_TEXT
        *
        results[
            "probability_roberta"
        ]
        +
        ALPHA_IMAGE
        *
        results[
            "probability_resnet"
        ]
    )


    results[
        "prediction_fusion"
    ] = (
        results[
            "probability_fusion"
        ]
        >= THRESHOLD
    ).astype(int)


    labels = (
        results[
            "label"
        ].to_numpy()
    )


    # ========================================================
    # Metrics
    # ========================================================

    systems = {
        "roberta": (
            results[
                "prediction_roberta"
            ].to_numpy(),

            results[
                "probability_roberta"
            ].to_numpy(),
        ),

        "resnet": (
            results[
                "prediction_resnet"
            ].to_numpy(),

            results[
                "probability_resnet"
            ].to_numpy(),
        ),

        "late_fusion": (
            results[
                "prediction_fusion"
            ].to_numpy(),

            results[
                "probability_fusion"
            ].to_numpy(),
        ),
    }


    metrics = {}


    print(
        "\n" + "=" * 70
    )

    print(
        "FINAL PERFORMANCE"
    )

    print("=" * 70)


    for name, (
        predictions,
        probabilities
    ) in systems.items():

        model_metrics = (
            calculate_metrics(
                labels,
                predictions,
                probabilities
            )
        )

        model_metrics[
            "ece"
        ] = (
            expected_calibration_error(
                labels,
                probabilities
            )
        )

        metrics[
            name
        ] = model_metrics


        print(
            "\n" + name.upper()
        )

        print(
            "-" * len(name)
        )


        for key in [
            "accuracy",
            "precision",
            "recall",
            "f1",
            "f1_macro",
            "roc_auc",
            "pr_auc",
            "brier_score",
            "log_loss",
            "ece",
        ]:

            print(
                f"{key:12s}: "
                f"{model_metrics[key]:.4f}"
            )


        print(
            "Confusion matrix:"
        )

        print(
            np.array(
                model_metrics[
                    "confusion_matrix"
                ]
            )
        )


    # ========================================================
    # Final paired significance:
    # late fusion vs RoBERTa
    # ========================================================

    roberta_pred = (
        systems[
            "roberta"
        ][0]
    )

    roberta_prob = (
        systems[
            "roberta"
        ][1]
    )

    fusion_pred = (
        systems[
            "late_fusion"
        ][0]
    )

    fusion_prob = (
        systems[
            "late_fusion"
        ][1]
    )


    roberta_correct = (
        roberta_pred
        == labels
    )

    fusion_correct = (
        fusion_pred
        == labels
    )


    roberta_only = int(
        np.sum(
            roberta_correct
            &
            ~fusion_correct
        )
    )

    fusion_only = int(
        np.sum(
            ~roberta_correct
            &
            fusion_correct
        )
    )


    discordant = (
        roberta_only
        +
        fusion_only
    )


    if discordant > 0:

        mcnemar_p = float(
            binomtest(
                min(
                    roberta_only,
                    fusion_only
                ),
                n=discordant,
                p=0.5,
                alternative="two-sided"
            ).pvalue
        )

    else:

        mcnemar_p = 1.0


    print(
        "\n" + "=" * 70
    )

    print(
        "FINAL FUSION VS ROBERTA "
        "PAIRED COMPARISON"
    )

    print("=" * 70)


    print(
        "\nRoBERTa correct / "
        "Fusion wrong:",
        roberta_only
    )

    print(
        "RoBERTa wrong / "
        "Fusion correct:",
        fusion_only
    )

    print(
        "Discordant:",
        discordant
    )

    print(
        f"McNemar exact p-value: "
        f"{mcnemar_p:.6f}"
    )


    observed_differences = {}


    print(
        "\nObserved differences "
        "(Fusion - RoBERTa):"
    )


    for metric in [
        "accuracy",
        "f1",
        "f1_macro",
        "roc_auc",
        "pr_auc",
    ]:

        difference = (
            metrics[
                "late_fusion"
            ][metric]
            -
            metrics[
                "roberta"
            ][metric]
        )

        observed_differences[
            metric
        ] = float(
            difference
        )

        print(
            f"{metric:12s}: "
            f"{difference:+.4f}"
        )


    print(
        f"\nRunning "
        f"{BOOTSTRAP_SAMPLES:,} "
        "paired bootstrap samples..."
    )


    bootstrap = paired_bootstrap(
        labels,
        roberta_pred,
        roberta_prob,
        fusion_pred,
        fusion_prob
    )


    print(
        "\n95% paired bootstrap "
        "confidence intervals:"
    )


    for metric in [
        "accuracy",
        "f1",
        "f1_macro",
        "roc_auc",
        "pr_auc",
    ]:

        lower = (
            bootstrap[
                metric
            ][
                "ci_95_lower"
            ]
        )

        upper = (
            bootstrap[
                metric
            ][
                "ci_95_upper"
            ]
        )

        observed = (
            observed_differences[
                metric
            ]
        )


        print(
            f"{metric:12s}: "
            f"{observed:+.4f} "
            f"[{lower:+.4f}, "
            f"{upper:+.4f}]"
        )


    # ========================================================
    # Save final outputs
    # ========================================================

    results.to_csv(
        OUTPUT_ROOT
        / "final_predictions.csv",
        index=False
    )


    final_output = {
        "holdout": {
            "samples":
                int(
                    len(results)
                ),

            "ordered_id_sha256":
                fingerprint,

            "label_counts": {
                str(key):
                    int(value)

                for key, value
                in dataframe[
                    "label"
                ]
                .value_counts()
                .sort_index()
                .items()
            },
        },

        "locked_specification": {
            "alpha_text":
                ALPHA_TEXT,

            "alpha_image":
                ALPHA_IMAGE,

            "threshold":
                THRESHOLD,

            "max_length":
                MAX_LENGTH,

            "image_size":
                224,
        },

        "metrics":
            metrics,

        "fusion_vs_roberta": {
            "roberta_correct_fusion_wrong":
                roberta_only,

            "roberta_wrong_fusion_correct":
                fusion_only,

            "discordant":
                discordant,

            "mcnemar_exact_p":
                mcnemar_p,

            "observed_differences":
                observed_differences,

            "bootstrap_samples":
                BOOTSTRAP_SAMPLES,

            "bootstrap_ci_95":
                bootstrap,
        },
    }


    with (
        OUTPUT_ROOT
        / "final_results.json"
    ).open(
        "w",
        encoding="utf-8"
    ) as f:

        json.dump(
            final_output,
            f,
            indent=2
        )


    print(
        "\n" + "=" * 70
    )

    print(
        "FINAL EVALUATION COMPLETE"
    )

    print("=" * 70)

    print(
        "\nResults saved to:",
        OUTPUT_ROOT
    )

    print(
        "\nThese are the locked final "
        "holdout results."
    )


# END REGISTERED SOURCE BLOCK


In [76]:
%%project_source multimodal-fake-news-detection/scripts/evaluate_final_holdout.py 4
if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


<a id="methodology"></a>
## 8. Later methodology notebook

The original explanatory Markdown and all eight code cells are reproduced below. They run as one separate notebook when explicitly requested, because later cells depend on earlier variables. The initial setup resolves the original-project and v2 folders relative to a repository root. Outputs and manifests are written under that working copy. Embedded original outputs are omitted; saved evidence is available separately below.

# Fakeddit multimodal methodology audit — v2

This notebook adds the methodological checks that were missing from the original project while preserving the original code, data, checkpoints, and results. It reads from the sibling `multimodal-fake-news-detection` folder and writes only to this `v2` folder.

The notebook covers:

1. binary-label semantics and internal consistency;
2. class-dependent image-selection bias;
3. a fairer validation-tuned and calibrated RoBERTa comparison;
4. source, domain, and time subgroup performance plus a source-only shortcut baseline;
5. perceptual-image duplicate screening;
6. source-disjoint and chronological manifests for stronger future retraining;
7. explainability coverage and reporting consistency checks.

The final holdout is used only for locked evaluation of predeclared controls. No original model or result is overwritten.

**Original methodology code cell 1**

In [77]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell1 0
from pathlib import Path
import json, hashlib, math, warnings
import numpy as np
import pandas as pd
import matplotlib.pyplot as plt
from PIL import Image
from scipy.fft import dctn
from scipy.stats import chi2_contingency
from sklearn.calibration import calibration_curve
from sklearn.linear_model import LogisticRegression
from sklearn.metrics import (
    accuracy_score, precision_score, recall_score, f1_score,
    roc_auc_score, average_precision_score, brier_score_loss,
    log_loss, confusion_matrix
)
from sklearn.model_selection import train_test_split

# Open the notebook from v2 or the submission repository root.
REPO_ROOT = Path.cwd().resolve()
if REPO_ROOT.name == "v2":
    REPO_ROOT = REPO_ROOT.parent
ORIGINAL_ROOT = REPO_ROOT / "multimodal-fake-news-detection"
V2_ROOT = REPO_ROOT / "v2"
OUTPUT_ROOT = V2_ROOT / "outputs"
MANIFEST_ROOT = V2_ROOT / "manifests"
RAW_ROOT = ORIGINAL_ROOT / "data" / "raw" / "fakeddit"
PROCESSED_ROOT = ORIGINAL_ROOT / "data" / "processed" / "fakeddit"
RESULTS_ROOT = ORIGINAL_ROOT / "results"
SEED = 2026

assert ORIGINAL_ROOT.exists(), ORIGINAL_ROOT
assert V2_ROOT != ORIGINAL_ROOT and ORIGINAL_ROOT not in V2_ROOT.parents
OUTPUT_ROOT.mkdir(parents=True, exist_ok=True)
MANIFEST_ROOT.mkdir(parents=True, exist_ok=True)

def save_json(name, obj):
    path = OUTPUT_ROOT / name
    path.write_text(json.dumps(obj, indent=2, default=str), encoding="utf-8")
    return path

def raw_path(split):
    name = {"train":"multimodal_train.tsv", "validation":"multimodal_validate.tsv", "test":"multimodal_test_public.tsv"}[split]
    return RAW_ROOT / "multimodal_only_samples" / name

def read_raw(split, columns=None):
    return pd.read_csv(raw_path(split), sep="\t", usecols=columns, low_memory=False)

def metrics(y, p, threshold=0.5):
    y = np.asarray(y, dtype=int); p = np.clip(np.asarray(p, dtype=float), 1e-7, 1-1e-7)
    pred = (p >= threshold).astype(int)
    return {
        "n": int(len(y)), "threshold": float(threshold),
        "accuracy": float(accuracy_score(y, pred)),
        "precision": float(precision_score(y, pred, zero_division=0)),
        "recall": float(recall_score(y, pred, zero_division=0)),
        "f1": float(f1_score(y, pred, zero_division=0)),
        "macro_f1": float(f1_score(y, pred, average="macro", zero_division=0)),
        "roc_auc": float(roc_auc_score(y, p)) if len(np.unique(y)) == 2 else np.nan,
        "pr_auc": float(average_precision_score(y, p)) if len(np.unique(y)) == 2 else np.nan,
        "brier": float(brier_score_loss(y, p)),
        "log_loss": float(log_loss(y, p, labels=[0,1])),
        "confusion_matrix": confusion_matrix(y, pred, labels=[0,1]).tolist(),
    }

print("Original (read-only):", ORIGINAL_ROOT)
print("v2 outputs:", V2_ROOT)
# END REGISTERED SOURCE BLOCK


## 1. Verify label semantics

Fakeddit's six-way label `0` is the true-content category; the other five categories are forms of false or misleading content. The binary encoding is therefore checked programmatically: binary class `1` must correspond exactly to six-way class `0`, and binary class `0` to six-way classes `1–5`.

**Original methodology code cell 3**

In [78]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell3 0
label_rows = []
label_tables = {}
for split in ["train", "validation", "test"]:
    d = read_raw(split, ["id", "2_way_label", "3_way_label", "6_way_label"])
    tab = pd.crosstab(d["2_way_label"], d["6_way_label"])
    label_tables[split] = tab
    consistent = ((d["2_way_label"] == 1) == (d["6_way_label"] == 0))
    label_rows.append({
        "split": split, "n": len(d), "consistent_n": int(consistent.sum()),
        "inconsistent_n": int((~consistent).sum()), "consistent_pct": float(100*consistent.mean())
    })
    display(tab)

label_audit = pd.DataFrame(label_rows)
label_audit.to_csv(OUTPUT_ROOT / "label_semantics_audit.csv", index=False)
assert label_audit["inconsistent_n"].sum() == 0
semantics = {
    "binary_class_1": "true/real content",
    "binary_class_0": "fake or misleading content (six-way classes 1-5)",
    "verification": label_rows,
    "limitation": "This verifies dataset encoding, not the factual correctness of every distant-supervision label."
}
save_json("label_semantics.json", semantics)
display(label_audit)
# END REGISTERED SOURCE BLOCK


## 2. Quantify selection bias caused by image availability

Equal sample IDs make comparisons between modalities fair within the retained subset. They do not make that subset representative. This section measures retention by label, year, domain, and subreddit and tests whether retention is independent of the binary label.

**Original methodology code cell 5**

In [79]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell5 0
status_parts = []
for split in ["train", "validation", "test"]:
    p = PROCESSED_ROOT / "development_clean" / f"{split}_with_image_status.parquet"
    s = pd.read_parquet(p)
    meta = read_raw(split, ["id", "subreddit", "domain", "created_utc", "2_way_label"])
    s["id"] = s["id"].astype(str); meta["id"] = meta["id"].astype(str)
    s = s.merge(meta, on="id", how="left", validate="one_to_one")
    s["retained"] = s["image_usable"].fillna(False).astype(bool)
    s["year"] = pd.to_datetime(s["created_utc"], unit="s", errors="coerce", utc=True).dt.year
    status_parts.append(s)
status = pd.concat(status_parts, ignore_index=True)

retention = (status.groupby(["split", "label"])["retained"]
             .agg(total="size", retained="sum", retention_rate="mean").reset_index())
retention["removed"] = retention["total"] - retention["retained"]
retention.to_csv(OUTPUT_ROOT / "selection_retention_by_label.csv", index=False)

contingency = pd.crosstab(status["label"], status["retained"])
chi2, p_value, _, _ = chi2_contingency(contingency)
n = contingency.to_numpy().sum()
cramers_v = math.sqrt(chi2 / n)
bias_summary = {
    "n": int(n), "chi_square": float(chi2), "p_value": float(p_value),
    "cramers_v": float(cramers_v),
    "interpretation": "Large dependence means complete-case filtering changes the target population. Macro-F1 does not remove this selection bias."
}
save_json("selection_bias_summary.json", bias_summary)

for group in ["subreddit", "domain", "year"]:
    g = (status.groupby(group, dropna=False)["retained"]
         .agg(total="size", retained="sum", retention_rate="mean").reset_index())
    g["removed"] = g["total"] - g["retained"]
    g.sort_values(["total", "retention_rate"], ascending=[False, True]).to_csv(
        OUTPUT_ROOT / f"selection_retention_by_{group}.csv", index=False)

display(retention)
print(bias_summary)

fig, ax = plt.subplots(figsize=(7,4))
for split, grp in retention.groupby("split"):
    ax.plot(grp["label"].astype(str), grp["retention_rate"], marker="o", label=split)
ax.set(xlabel="Binary label (0=fake/misleading, 1=true)", ylabel="Image retention rate", ylim=(0,1),
       title="Image filtering is strongly class-dependent")
ax.legend(); fig.tight_layout()
fig.savefig(OUTPUT_ROOT / "selection_retention_by_label.png", dpi=180)
plt.show()
# END REGISTERED SOURCE BLOCK


## 3. Fair text-only threshold and calibration controls

The original fusion weight was selected on validation macro-F1 while RoBERTa used the default 0.5 threshold. This section gives RoBERTa the same opportunity to tune its decision threshold. It also fits Platt calibration on one stratified half of validation and selects its threshold on the other half, then evaluates each predeclared variant once on the frozen holdout.

**Original methodology code cell 7**

In [80]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell7 0
val = pd.read_csv(RESULTS_ROOT / "metrics" / "baseline_probabilities" / "roberta_validation.csv")
final = pd.read_csv(RESULTS_ROOT / "metrics" / "final_evaluation" / "final_predictions.csv")
val = val.rename(columns={"probability_class_1":"p_text"})

threshold_grid = np.linspace(0.05, 0.95, 181)
threshold_scores = pd.DataFrame({
    "threshold": threshold_grid,
    "validation_macro_f1": [metrics(val.label, val.p_text, t)["macro_f1"] for t in threshold_grid]
})
best_t = float(threshold_scores.sort_values(["validation_macro_f1", "threshold"], ascending=[False, True]).iloc[0].threshold)
threshold_scores.to_csv(OUTPUT_ROOT / "roberta_validation_threshold_search.csv", index=False)

idx_cal, idx_tune = train_test_split(np.arange(len(val)), test_size=0.5, random_state=SEED, stratify=val.label)
def logit(p):
    p = np.clip(np.asarray(p, float), 1e-6, 1-1e-6)
    return np.log(p/(1-p)).reshape(-1,1)
platt = LogisticRegression(C=1e6, solver="lbfgs", random_state=SEED)
platt.fit(logit(val.p_text.iloc[idx_cal]), val.label.iloc[idx_cal])
p_tune = platt.predict_proba(logit(val.p_text.iloc[idx_tune]))[:,1]
platt_grid = pd.DataFrame({
    "threshold": threshold_grid,
    "tuning_half_macro_f1": [metrics(val.label.iloc[idx_tune], p_tune, t)["macro_f1"] for t in threshold_grid]
})
platt_t = float(platt_grid.sort_values(["tuning_half_macro_f1", "threshold"], ascending=[False, True]).iloc[0].threshold)
platt_grid.to_csv(OUTPUT_ROOT / "roberta_platt_threshold_search.csv", index=False)
p_final_platt = platt.predict_proba(logit(final.probability_roberta))[:,1]

control_results = {
    "roberta_default_0.5": metrics(final.label, final.probability_roberta, 0.5),
    "roberta_validation_tuned_threshold": metrics(final.label, final.probability_roberta, best_t),
    "roberta_platt_default_0.5": metrics(final.label, p_final_platt, 0.5),
    "roberta_platt_tuned_threshold": metrics(final.label, p_final_platt, platt_t),
    "locked_late_fusion": metrics(final.label, final.probability_fusion, 0.5),
}
control_table = pd.DataFrame(control_results).T.reset_index(names="model")
control_table.to_csv(OUTPUT_ROOT / "fair_text_baseline_comparison.csv", index=False)
save_json("fair_text_baseline_comparison.json", {
    "validation_selected_text_threshold": best_t,
    "platt_calibration_fit_n": int(len(idx_cal)), "platt_threshold_tuning_n": int(len(idx_tune)),
    "platt_selected_threshold": platt_t, "final_results": control_results
})
display(control_table[["model","accuracy","macro_f1","roc_auc","pr_auc","brier","log_loss","threshold"]])
# END REGISTERED SOURCE BLOCK


## 4. Source, domain, and time diagnostics

These are subgroup diagnostics, not a source-disjoint test: the trained models may have seen the same source categories during training. A source-only baseline is also fitted from original training labels. If it performs well, source identity alone carries target information and remains a plausible shortcut even though metadata was withheld from the neural networks.

**Original methodology code cell 9**

In [81]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell9 0
test_meta = read_raw("test", ["id","subreddit","domain","created_utc","2_way_label"])
test_meta["id"] = test_meta["id"].astype(str); final["id"] = final["id"].astype(str)
enriched = final.merge(test_meta, on="id", how="left", validate="one_to_one")
enriched["year"] = pd.to_datetime(enriched.created_utc, unit="s", errors="coerce", utc=True).dt.year

def subgroup_table(group, min_n=30):
    rows=[]
    for key, g in enriched.groupby(group, dropna=False):
        if len(g) < min_n or g.label.nunique() < 2: continue
        tm=metrics(g.label, g.probability_roberta); fm=metrics(g.label, g.probability_fusion)
        rows.append({group:key, "n":len(g), "class_1_rate":g.label.mean(),
                     "roberta_macro_f1":tm["macro_f1"], "fusion_macro_f1":fm["macro_f1"],
                     "fusion_delta_macro_f1":fm["macro_f1"]-tm["macro_f1"],
                     "roberta_accuracy":tm["accuracy"], "fusion_accuracy":fm["accuracy"]})
    columns=[group,"n","class_1_rate","roberta_macro_f1","fusion_macro_f1",
             "fusion_delta_macro_f1","roberta_accuracy","fusion_accuracy"]
    return pd.DataFrame(rows, columns=columns).sort_values("n", ascending=False)

for group in ["subreddit","domain","year"]:
    table=subgroup_table(group)
    table.to_csv(OUTPUT_ROOT / f"final_performance_by_{group}.csv", index=False)
    display(table.head(15))

train_source = read_raw("train", ["subreddit","2_way_label"])
global_rate = float(train_source["2_way_label"].mean())
rates = train_source.groupby("subreddit")["2_way_label"].agg(["mean","size"])
smooth = (rates["mean"]*rates["size"] + global_rate*50)/(rates["size"]+50)
source_prob = enriched["subreddit"].map(smooth).fillna(global_rate).to_numpy()
source_only = metrics(enriched.label, source_prob, 0.5)

source_label_tab = pd.crosstab(train_source.subreddit, train_source["2_way_label"])
chi2, p, _, _ = chi2_contingency(source_label_tab)
v = math.sqrt(chi2/(source_label_tab.to_numpy().sum()*min(source_label_tab.shape[0]-1, source_label_tab.shape[1]-1)))
source_summary={"source_only_final_holdout":source_only,"training_source_label_cramers_v":float(v),"chi_square_p":float(p)}
save_json("source_shortcut_audit.json", source_summary)
print(source_summary)
# END REGISTERED SOURCE BLOCK


## 5. Perceptual duplicate screening

Exact hashes miss resized or recompressed copies. A 64-bit perceptual hash is computed for every usable development image and final image. A BK-tree searches for cross-set pairs within Hamming distance 6. These pairs are candidates for manual review; perceptual similarity alone is not proof of duplication.

**Original methodology code cell 11**

In [82]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell11 0
def resolve_original(path_value):
    p=Path(str(path_value)); return p if p.is_absolute() else ORIGINAL_ROOT/p

def phash64(path):
    with Image.open(path) as im:
        a=np.asarray(im.convert("L").resize((32,32), Image.Resampling.LANCZOS), dtype=float)
    low=dctn(a, type=2, norm="ortho")[:8,:8]
    med=np.median(low.ravel()[1:])
    bits=(low>med).ravel()
    value=0
    for bit in bits: value=(value<<1)|int(bit)
    return value

cache_path=OUTPUT_ROOT/"perceptual_hashes.csv"
if cache_path.exists():
    hashes=pd.read_csv(cache_path, dtype={"id":str,"phash_hex":str})
else:
    image_rows=[]
    for split in ["train","validation","test"]:
        d=pd.read_parquet(PROCESSED_ROOT/"development_clean"/f"{split}.parquet")
        image_rows.extend(("development",str(r.id),resolve_original(r.image_path)) for r in d.itertuples())
    hold=pd.read_parquet(PROCESSED_ROOT/"final_holdout"/"final_5000.parquet")
    image_rows.extend(("final",str(r.id),resolve_original(r.image_path)) for r in hold.itertuples())
    out=[]
    for i,(partition,sid,path) in enumerate(image_rows,1):
        try: out.append({"partition":partition,"id":sid,"path":str(path),"phash_hex":f"{phash64(path):016x}","error":""})
        except Exception as e: out.append({"partition":partition,"id":sid,"path":str(path),"phash_hex":"","error":type(e).__name__})
        if i%2500==0: print(f"Hashed {i:,}/{len(image_rows):,}")
    hashes=pd.DataFrame(out); hashes.to_csv(cache_path,index=False)

class BKNode:
    def __init__(self,key,payload): self.key,self.payload,self.children=key,[payload],{}
    def add(self,key,payload):
        node=self
        while True:
            dist=(node.key^key).bit_count()
            if dist==0: node.payload.append(payload); return
            if dist not in node.children: node.children[dist]=BKNode(key,payload); return
            node=node.children[dist]
    def search(self,key,radius):
        found=[]; stack=[self]
        while stack:
            node=stack.pop(); dist=(node.key^key).bit_count()
            if dist<=radius: found.extend((p,dist) for p in node.payload)
            stack.extend(child for edge,child in node.children.items() if dist-radius<=edge<=dist+radius)
        return found

dev=hashes[(hashes.partition=="development") & hashes.phash_hex.ne("")]
fin=hashes[(hashes.partition=="final") & hashes.phash_hex.ne("")]
tree=None
for r in dev.itertuples():
    key=int(r.phash_hex,16)
    if tree is None: tree=BKNode(key,(r.id,r.path,r.phash_hex))
    else: tree.add(key,(r.id,r.path,r.phash_hex))
pairs=[]
for r in fin.itertuples():
    for (dev_id,dev_path,dev_hash),distance in tree.search(int(r.phash_hex,16),6):
        pairs.append({"final_id":r.id,"development_id":dev_id,"hamming_distance":distance,
                      "final_path":r.path,"development_path":dev_path,"final_phash":r.phash_hex,"development_phash":dev_hash})
near=pd.DataFrame(pairs).sort_values(["hamming_distance","final_id"]) if pairs else pd.DataFrame(columns=["final_id","development_id","hamming_distance"])
near.to_csv(OUTPUT_ROOT/"perceptual_near_duplicate_candidates.csv",index=False)
print(f"Usable hashes: development={len(dev):,}; final={len(fin):,}")
print(f"Cross-set candidate pairs at Hamming distance <=6: {len(near):,}")
display(near.head(20))
# END REGISTERED SOURCE BLOCK


## 6. Stronger split manifests for future retraining

The current checkpoints cannot be converted into source-disjoint or chronological experiments after training. This section creates reproducible manifests for those experiments without running expensive model training. Each manifest uses only the existing cleaned multimodal development examples.

**Original methodology code cell 13**

In [83]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell13 0
clean_parts=[]
for split in ["train","validation","test"]:
    d=pd.read_parquet(PROCESSED_ROOT/"development_clean"/f"{split}.parquet")
    meta=read_raw(split,["id","subreddit","domain","created_utc","2_way_label"])
    d["id"]=d.id.astype(str); meta["id"]=meta.id.astype(str)
    clean_parts.append(d.merge(meta,on="id",how="left",validate="one_to_one"))
clean=pd.concat(clean_parts,ignore_index=True).drop_duplicates("id")
clean["created_datetime"]=pd.to_datetime(clean.created_utc,unit="s",errors="coerce",utc=True)

# Source-disjoint: Fakeddit subreddits are label-pure. Allocate whole subreddits
# separately inside each label so every split contains both classes.
purity=clean.groupby("subreddit")["label"].nunique()
assert purity.max()==1, "Expected subreddit-level distant-supervision labels."
source_labels=clean.groupby("subreddit")["label"].first()
counts=clean.groupby("subreddit").size()
assignment={}
for label in sorted(clean.label.unique()):
    label_counts=counts[source_labels==label].sort_values(ascending=False)
    label_total=int(label_counts.sum())
    targets={"train":.70*label_total,"validation":.15*label_total,"test":.15*label_total}
    totals={k:0 for k in targets}
    for source,count in label_counts.items():
        split=min(targets,key=lambda k: totals[k]/targets[k])
        assignment[source]=split; totals[split]+=int(count)
source_manifest=clean[["id","label","text","image_path","subreddit","domain","created_utc"]].copy()
source_manifest["v2_split"]=source_manifest.subreddit.map(assignment)
assert source_manifest.groupby("subreddit").v2_split.nunique().max()==1
assert source_manifest.groupby("v2_split").label.nunique().min()==2
source_manifest.to_parquet(MANIFEST_ROOT/"source_disjoint.parquet",index=False)

chronological=clean.sort_values(["created_datetime","id"]).copy()
chronological["v2_split"]="train"
chronological.iloc[int(.70*len(chronological)):int(.85*len(chronological)), chronological.columns.get_loc("v2_split")]="validation"
chronological.iloc[int(.85*len(chronological)):, chronological.columns.get_loc("v2_split")]="test"
chronological[["id","label","text","image_path","subreddit","domain","created_utc","v2_split"]].to_parquet(
    MANIFEST_ROOT/"chronological.parquet",index=False)

split_summary=pd.concat([
    source_manifest.groupby("v2_split").agg(n=("id","size"),class_1_rate=("label","mean")).assign(manifest="source_disjoint"),
    chronological.groupby("v2_split").agg(n=("id","size"),class_1_rate=("label","mean")).assign(manifest="chronological")
]).reset_index()
split_summary.to_csv(OUTPUT_ROOT/"v2_manifest_summary.csv",index=False)
display(split_summary)
# END REGISTERED SOURCE BLOCK


## 7. Explainability coverage and reporting checks

This verifies whether the stored artifacts match the method description and writes a machine-readable correction list for the dissertation draft.

**Original methodology code cell 15**

In [84]:
%%project_source v2/methodology_gap_analysis_v2.ipynb::cell15 0
cases32=pd.read_csv(RESULTS_ROOT/"case_studies"/"all_32_multimodal_cases.csv")
cases8=pd.read_csv(RESULTS_ROOT/"case_studies"/"selected_8_case_studies.csv")
shap_summary=pd.read_csv(RESULTS_ROOT/"shap"/"shap_case_summary.csv")
grad_summary=pd.read_csv(RESULTS_ROOT/"gradcam"/"gradcam_case_summary.csv")
coverage={
    "all_multimodal_cases":int(len(cases32)), "selected_paired_cases":int(len(cases8)),
    "shap_cases":int(len(shap_summary)), "gradcam_cases":int(len(grad_summary)),
    "case_columns":list(cases32.columns),
}
if "label" in cases32.columns: coverage["all_32_label_counts"]={str(k):int(v) for k,v in cases32.label.value_counts().items()}
save_json("explainability_coverage.json",coverage)

raw_test_n=len(read_raw("test",["id"]))
robustness=json.loads((RESULTS_ROOT/"metrics"/"missing_modality_robustness"/"results.json").read_text())
changes={r["scenario"]:r["macro_f1_change_vs_full"] for r in robustness["results"]}
checks=pd.DataFrame([
    {"item":"public test size","observed":raw_test_n,"expected":59319,"status":"PASS" if raw_test_n==59319 else "FAIL","draft_action":"Use 59,319 consistently."},
    {"item":"missing text change sign","observed":changes.get("missing_text_image_fallback"),"expected":"negative","status":"PASS" if changes.get("missing_text_image_fallback",1)<0 else "FAIL","draft_action":"Report -0.0906, not +0.0906."},
    {"item":"32-case table exists","observed":len(cases32),"expected":32,"status":"PASS" if len(cases32)==32 else "FAIL","draft_action":"Describe the full 32-case analysis and distinguish it from the four illustrated cases."},
    {"item":"paired SHAP and Grad-CAM coverage","observed":f"SHAP={len(shap_summary)}, Grad-CAM={len(grad_summary)}","expected":">=32 each","status":"PASS" if min(len(shap_summary),len(grad_summary))>=32 else "FAIL","draft_action":"Reconcile claimed and generated explanation counts."},
])
checks.to_csv(OUTPUT_ROOT/"reporting_consistency_checks.csv",index=False)
display(checks)
print(coverage)
# END REGISTERED SOURCE BLOCK


## Interpretation boundaries

The strongest supported conclusion remains specific: on the selected cleaned Fakeddit sample and locked checkpoints, late probability fusion improves over the original RoBERTa decision rule. The added controls show whether that advantage remains after fair threshold tuning and how strongly source and selection effects constrain generalisation.

The source-disjoint and chronological manifests must be used to retrain all models from scratch before making claims about transfer to unseen sources or later periods. Full training-seed uncertainty likewise requires several independent end-to-end training runs; it cannot be recovered from one checkpoint. This notebook deliberately does not fabricate those results.

<a id="source"></a>
## 9. Source-disjoint retraining

This runner implements `audit â†’ smoke â†’ train-roberta â†’ train-resnet â†’ lock â†’ test`. Both encoders are retrained on the new training partition. The validation partition determines the coefficient, even when its choice later performs poorly on test. The submission version replaces hard-coded original paths with repository-relative paths and an optional `FAKEDDIT_PROJECT_ROOT`; the earlier local version is preserved in the appendix.

### 9.1 Run source disjoint

Audit the source-disjoint manifests, smoke-test inputs, retrain both encoders, lock fusion on validation and evaluate the separate test partition.

**Source:** `v2/experiments/source_disjoint/run_source_disjoint.py`  
**Imported modules:** `PIL`, `__future__`, `argparse`, `datetime`, `hashlib`, `json`, `matplotlib`, `numpy`, `os`, `pandas`, `pathlib`, `platform`, `random`, `scipy`, `shutil`, `sklearn`, `sys`, `torch`, `torchvision`, `transformers`  
**Top-level components:** `paths`, `make_dirs`, `dump_json`, `set_seed`, `resolve_image_path`, `load_manifest`, `split_df`, `metrics_for`, `TextDataset`, `ImageDataset`, `image_transform`, `worker_seed`, `text_evaluate`, `image_evaluate`, `prediction_frame`, `stage_audit`, `create_resnet`, `stage_smoke`, `train_roberta`, `train_resnet`, `stage_lock`, `ece`, `calibration_for`, `bootstrap`, `reliability_plot`, `markdown_table`, `stage_test`, `main`

The following cells contain the complete source; Run All registers it for inspection/export.

In [85]:
%%project_source v2/experiments/source_disjoint/run_source_disjoint.py 0
"""Isolated source-disjoint retraining and evaluation for the Fakeddit study.

The command is deliberately split into stages so the test partition is not used
until both validation checkpoints and the late-fusion coefficient are locked.
"""

from __future__ import annotations

import argparse
import hashlib
import json
import os
import platform
import random
import shutil
import sys
from datetime import datetime, timezone
from pathlib import Path

import matplotlib.pyplot as plt
import numpy as np
import pandas as pd
import scipy
import sklearn
import torch
import torch.nn as nn
import torchvision
import transformers
from PIL import Image
from scipy.stats import binomtest
from sklearn.linear_model import LogisticRegression
from sklearn.metrics import (
    accuracy_score,
    average_precision_score,
    brier_score_loss,
    confusion_matrix,
    f1_score,
    log_loss,
    precision_score,
    recall_score,
    roc_auc_score,
)
from torch.optim import AdamW
from torch.utils.data import DataLoader, Dataset
from torchvision import transforms
from torchvision.models import ResNet50_Weights, resnet50
from transformers import (
    AutoModelForSequenceClassification,
    AutoTokenizer,
    get_linear_schedule_with_warmup,
)


SEED = 42
MODEL_NAME = "roberta-base"
MAX_LENGTH = 64
THRESHOLD = 0.50
N_BINS = 10
N_BOOTSTRAPS = 5000
PLACEHOLDER_SHA256 = "faa24ec881e6040655c187a681d6dc496eb8aa41e1bd0652a180b3a40b457187"
REPOSITORY_ROOT = Path(__file__).resolve().parents[3]
PROJECT_ROOT = Path(os.environ.get("FAKEDDIT_PROJECT_ROOT", str(REPOSITORY_ROOT / "multimodal-fake-news-detection")))
SOURCE_MANIFEST = REPOSITORY_ROOT / "v2" / "manifests" / "source_disjoint.parquet"
DEFAULT_EXPERIMENT_ROOT = Path(__file__).resolve().parent


def paths(root: Path) -> dict[str, Path]:
    return {
        "root": root,
        "manifests": root / "manifests",
        "checkpoints": root / "checkpoints",
        "roberta_checkpoint": root / "checkpoints" / "roberta",
        "resnet_checkpoint": root / "checkpoints" / "resnet50",
        "predictions": root / "predictions",
        "metrics": root / "metrics",
        "logs": root / "logs",
        "figures": root / "figures",
        "bootstrap": root / "bootstrap",
        "calibration": root / "calibration",
        "reports": root / "reports",
        "manifest": root / "manifests" / "source_disjoint.parquet",
        "config": root / "experiment_config.json",
        "audit": root / "manifests" / "manifest_audit.json",
        "lock": root / "metrics" / "validation_lock.json",
    }


def make_dirs(root: Path) -> None:
    for key, value in paths(root).items():
        if key not in {"manifest", "config", "audit", "lock"}:
            value.mkdir(parents=True, exist_ok=True)


def dump_json(path: Path, value: dict) -> None:
    path.parent.mkdir(parents=True, exist_ok=True)
    path.write_text(json.dumps(value, indent=2, allow_nan=False), encoding="utf-8")


def set_seed(seed: int = SEED) -> None:
    os.environ["PYTHONHASHSEED"] = str(seed)
    random.seed(seed)
    np.random.seed(seed)
    torch.manual_seed(seed)
    if torch.cuda.is_available():
        torch.cuda.manual_seed_all(seed)
    torch.backends.cudnn.deterministic = True
    torch.backends.cudnn.benchmark = False


def resolve_image_path(value: str) -> Path:
    # Archived manifests retain the original workstation's absolute image paths.
    normalised = str(value).replace("\\", "/")
    marker = "/multimodal-fake-news-detection/"
    if marker in normalised:
        return PROJECT_ROOT / normalised.split(marker, 1)[1]
    path = Path(normalised)
    return path if path.is_absolute() else PROJECT_ROOT / path


def load_manifest(root: Path) -> pd.DataFrame:
    path = paths(root)["manifest"]
    if not path.exists():
        raise FileNotFoundError(f"Run the audit stage first: {path}")
    df = pd.read_parquet(path)
    required = {"id", "label", "text", "image_path", "subreddit", "v2_split"}
    missing = required.difference(df.columns)
    if missing:
        raise ValueError(f"Manifest lacks columns: {sorted(missing)}")
    df = df.copy()
    df["id"] = df["id"].astype(str)
    df["label"] = df["label"].astype(int)
    df["resolved_image_path"] = df["image_path"].map(lambda x: str(resolve_image_path(x)))
    return df


def split_df(df: pd.DataFrame, split: str) -> pd.DataFrame:
    result = df.loc[df["v2_split"].eq(split)].copy().reset_index(drop=True)
    if result.empty:
        raise ValueError(f"Empty split: {split}")
    return result


def metrics_for(labels, predictions, probabilities) -> dict:
    labels = np.asarray(labels, dtype=int)
    predictions = np.asarray(predictions, dtype=int)
    probabilities = np.asarray(probabilities, dtype=float)
    result = {
        "accuracy": float(accuracy_score(labels, predictions)),
        "precision": float(precision_score(labels, predictions, zero_division=0)),
        "recall": float(recall_score(labels, predictions, zero_division=0)),
        "f1": float(f1_score(labels, predictions, zero_division=0)),
        "macro_f1": float(f1_score(labels, predictions, average="macro", zero_division=0)),
        "recall_class_0": float(recall_score(labels, predictions, labels=[0], average=None, zero_division=0)[0]),
        "recall_class_1": float(recall_score(labels, predictions, labels=[1], average=None, zero_division=0)[0]),
        "roc_auc": float(roc_auc_score(labels, probabilities)) if np.unique(labels).size == 2 else None,
        "pr_auc": float(average_precision_score(labels, probabilities)) if np.unique(labels).size == 2 else None,
        "confusion_matrix": confusion_matrix(labels, predictions, labels=[0, 1]).tolist(),
    }
    return result


# END REGISTERED SOURCE BLOCK


In [86]:
%%project_source v2/experiments/source_disjoint/run_source_disjoint.py 1
class TextDataset(Dataset):
    def __init__(self, dataframe: pd.DataFrame, tokenizer):
        self.ids = dataframe["id"].astype(str).tolist()
        self.labels = torch.tensor(dataframe["label"].to_numpy(dtype=int), dtype=torch.long)
        self.encodings = tokenizer(
            dataframe["text"].fillna("").astype(str).tolist(),
            padding="max_length",
            truncation=True,
            max_length=MAX_LENGTH,
            return_tensors="pt",
        )

    def __len__(self):
        return len(self.labels)

    def __getitem__(self, index):
        item = {key: value[index] for key, value in self.encodings.items()}
        item["labels"] = self.labels[index]
        item["sample_index"] = torch.tensor(index, dtype=torch.long)
        return item


class ImageDataset(Dataset):
    def __init__(self, dataframe: pd.DataFrame, transform):
        self.df = dataframe.reset_index(drop=True)
        self.transform = transform

    def __len__(self):
        return len(self.df)

    def __getitem__(self, index):
        row = self.df.iloc[index]
        with Image.open(row["resolved_image_path"]) as image:
            tensor = self.transform(image.convert("RGB"))
        return {
            "image": tensor,
            "label": torch.tensor(int(row["label"]), dtype=torch.long),
            "sample_index": torch.tensor(index, dtype=torch.long),
        }


def image_transform():
    return transforms.Compose([
        transforms.Resize((224, 224)),
        transforms.ToTensor(),
        transforms.Normalize(mean=[0.485, 0.456, 0.406], std=[0.229, 0.224, 0.225]),
    ])


def worker_seed(worker_id: int) -> None:
    worker_seed_value = SEED + worker_id
    np.random.seed(worker_seed_value)
    random.seed(worker_seed_value)


def text_evaluate(model, loader, device):
    model.eval()
    labels, predictions, probabilities, indices = [], [], [], []
    total_loss = 0.0
    with torch.no_grad():
        for batch in loader:
            index = batch.pop("sample_index")
            cpu_labels = batch["labels"].numpy()
            batch = {key: value.to(device, non_blocking=True) for key, value in batch.items()}
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                output = model(**batch)
            probability = torch.softmax(output.logits, dim=1)[:, 1]
            prediction = (probability >= THRESHOLD).long()
            total_loss += float(output.loss.item())
            indices.extend(index.numpy().tolist())
            labels.extend(cpu_labels.tolist())
            predictions.extend(prediction.cpu().numpy().tolist())
            probabilities.extend(probability.cpu().float().numpy().tolist())
    result = metrics_for(labels, predictions, probabilities)
    result["loss"] = total_loss / len(loader)
    return result, np.asarray(indices), np.asarray(labels), np.asarray(predictions), np.asarray(probabilities)


def image_evaluate(model, loader, device):
    model.eval()
    labels, predictions, probabilities, indices = [], [], [], []
    total_loss = 0.0
    criterion = nn.CrossEntropyLoss()
    with torch.no_grad():
        for batch in loader:
            image = batch["image"].to(device, non_blocking=True)
            label = batch["label"].to(device, non_blocking=True)
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                logits = model(image)
                loss = criterion(logits, label)
            probability = torch.softmax(logits, dim=1)[:, 1]
            prediction = (probability >= THRESHOLD).long()
            total_loss += float(loss.item())
            indices.extend(batch["sample_index"].numpy().tolist())
            labels.extend(label.cpu().numpy().tolist())
            predictions.extend(prediction.cpu().numpy().tolist())
            probabilities.extend(probability.cpu().float().numpy().tolist())
    result = metrics_for(labels, predictions, probabilities)
    result["loss"] = total_loss / len(loader)
    return result, np.asarray(indices), np.asarray(labels), np.asarray(predictions), np.asarray(probabilities)


def prediction_frame(dataframe, indices, labels, predictions, probabilities, prefix: str) -> pd.DataFrame:
    indexed = dataframe.iloc[indices].reset_index(drop=True)
    if not np.array_equal(indexed["label"].to_numpy(dtype=int), labels):
        raise ValueError(f"Label alignment failed for {prefix}")
    return pd.DataFrame({
        "sample_id": indexed["id"].astype(str),
        "true_label": labels,
        f"{prefix}_probability_class1": probabilities,
        f"{prefix}_prediction": predictions,
    })


def stage_audit(root: Path) -> None:
    make_dirs(root)
    p = paths(root)
    if not SOURCE_MANIFEST.exists():
        raise FileNotFoundError(SOURCE_MANIFEST)
    if p["manifest"].exists():
        if hashlib.sha256(p["manifest"].read_bytes()).hexdigest() != hashlib.sha256(SOURCE_MANIFEST.read_bytes()).hexdigest():
            raise FileExistsError(f"An unrelated manifest already exists at {p['manifest']}")
    else:
        shutil.copy2(SOURCE_MANIFEST, p["manifest"])

    df = pd.read_parquet(p["manifest"])
    required = ["id", "label", "text", "image_path", "subreddit", "domain", "created_utc", "v2_split"]
    if list(df.columns) != required:
        raise ValueError(f"Unexpected schema: {df.columns.tolist()}")
    if df["id"].astype(str).duplicated().any():
        raise ValueError("Duplicate sample IDs")
    if set(df["v2_split"]) != {"train", "validation", "test"}:
        raise ValueError("Unexpected split labels")
    if set(df["label"].astype(int)) != {0, 1}:
        raise ValueError("Unexpected class labels")

    source_sets = {name: set(group["subreddit"].astype(str)) for name, group in df.groupby("v2_split")}
    overlap = {}
    names = sorted(source_sets)
    for i, left in enumerate(names):
        for right in names[i + 1:]:
            overlap[f"{left}__{right}"] = sorted(source_sets[left] & source_sets[right])
    if any(overlap.values()):
        raise ValueError(f"Source overlap found: {overlap}")

    records, unreadable, placeholders = [], [], []
    for row in df.itertuples(index=False):
        image_path = resolve_image_path(row.image_path)
        exists = image_path.is_file()
        readable = False
        digest = None
        error = None
        if exists:
            try:
                with Image.open(image_path) as image:
                    image.verify()
                readable = True
                digest = hashlib.sha256(image_path.read_bytes()).hexdigest()
            except Exception as exc:  # recorded in audit output
                error = repr(exc)
        if not readable:
            unreadable.append({"id": str(row.id), "path": str(image_path), "error": error or "missing"})
        if digest == PLACEHOLDER_SHA256:
            placeholders.append(str(row.id))
        records.append({"v2_split": row.v2_split, "label": int(row.label), "readable": readable})
    checks = pd.DataFrame(records)
    split_rows = []
    for split in ["train", "validation", "test"]:
        part = df[df["v2_split"].eq(split)]
        verified = checks[checks["v2_split"].eq(split)]
        split_rows.append({
            "split": split,
            "manifest_samples": int(len(part)),
            "retained_samples": int(verified["readable"].sum()),
            "removed_samples": int((~verified["readable"]).sum()),
            "removed_class_0": 0,
            "removed_class_1": 0,
            "class_0": int(part["label"].eq(0).sum()),
            "class_1": int(part["label"].eq(1).sum()),
            "class_1_rate": float(part["label"].mean()),
            "sources": int(part["subreddit"].nunique()),
        })
    if unreadable or placeholders:
        raise ValueError(f"Manifest contains {len(unreadable)} unreadable and {len(placeholders)} placeholder images")
    pd.DataFrame(split_rows).to_csv(p["manifests"] / "split_counts.csv", index=False)

    manifest_sha = hashlib.sha256(p["manifest"].read_bytes()).hexdigest()
    audit = {
        "source_manifest": str(SOURCE_MANIFEST),
        "isolated_manifest": str(p["manifest"]),
        "sha256": manifest_sha,
        "schema": {column: str(dtype) for column, dtype in df.dtypes.items()},
        "rows": int(len(df)),
        "duplicate_ids": 0,
        "blank_text": int(df["text"].fillna("").astype(str).str.strip().eq("").sum()),
        "source_overlap": overlap,
        "unreadable_images": unreadable,
        "known_placeholder_images": placeholders,
        "splits": split_rows,
        "positive_class": "1 (true)",
        "negative_class": "0 (fake or misleading)",
        "note": "The manifest was constructed from the existing cleaned multimodal pool, so its manifest and retained counts are equal.",
    }
    dump_json(p["audit"], audit)
    config = {
        "experiment": "source_disjoint",
        "created_utc": datetime.now(timezone.utc).isoformat(),
        "seed": SEED,
        "project_root": str(PROJECT_ROOT),
        "source_manifest": str(SOURCE_MANIFEST),
        "isolated_manifest": str(p["manifest"]),
        "manifest_sha256": manifest_sha,
        "split_counts": {row["split"]: row["retained_samples"] for row in split_rows},
        "positive_class": 1,
        "classification_threshold": THRESHOLD,
        "roberta": {"base_model": MODEL_NAME, "pretrained_base_weights": True, "max_length": MAX_LENGTH, "batch_size": 16, "optimizer": "AdamW", "learning_rate": 2e-5, "weight_decay": 0.01, "gradient_clipping": 1.0, "warmup_fraction": 0.10, "max_epochs": 3, "selection_metric": "validation_macro_f1", "checkpoint": str(p["roberta_checkpoint"])},
        "resnet50": {"base_model": "resnet50", "weights": "IMAGENET1K_V2", "fine_tune": "full network", "input_size": [224, 224], "batch_size": 32, "optimizer": "AdamW", "learning_rate": 1e-4, "weight_decay": 0.01, "max_epochs": 3, "selection_metric": "validation_macro_f1", "checkpoint": str(p["resnet_checkpoint"] / "best_model.pt")},
        "fusion": {"formula": "alpha * p_text + (1 - alpha) * p_image", "alpha_search": [round(x, 2) for x in np.arange(0, 1.0001, 0.05)], "selection_metric": "validation_macro_f1", "tie_break": "closest to 0.50, then lower alpha", "selected_alpha": None},
        "calibration": {"ece_bins": N_BINS, "convention": "confidence bins from 0.5 to 1.0"},
        "bootstrap": {"iterations": N_BOOTSTRAPS, "seed": SEED, "paired": True},
        "packages": {"python": platform.python_version(), "torch": torch.__version__, "torchvision": torchvision.__version__, "transformers": transformers.__version__, "pandas": pd.__version__, "numpy": np.__version__, "scikit_learn": sklearn.__version__, "scipy": scipy.__version__},
        "hardware": {"cuda_available": torch.cuda.is_available(), "cuda_version": torch.version.cuda, "gpu": torch.cuda.get_device_name(0) if torch.cuda.is_available() else None},
    }
    dump_json(p["config"], config)
    print(pd.DataFrame(split_rows).to_string(index=False))
    print(f"Audit saved: {p['audit']}")


# END REGISTERED SOURCE BLOCK


In [87]:
%%project_source v2/experiments/source_disjoint/run_source_disjoint.py 2
def create_resnet() -> nn.Module:
    model = resnet50(weights=ResNet50_Weights.IMAGENET1K_V2)
    model.fc = nn.Linear(model.fc.in_features, 2)
    return model


def stage_smoke(root: Path) -> None:
    set_seed()
    df = load_manifest(root)
    train = split_df(df, "train").sample(n=32, random_state=SEED).reset_index(drop=True)
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    tokenizer = AutoTokenizer.from_pretrained(MODEL_NAME)
    text_loader = DataLoader(TextDataset(train, tokenizer), batch_size=8, shuffle=False)
    text_model = AutoModelForSequenceClassification.from_pretrained(MODEL_NAME, num_labels=2).to(device)
    text_batch = next(iter(text_loader))
    text_indices = text_batch.pop("sample_index")
    with torch.no_grad(), torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
        text_out = text_model(**{key: value.to(device) for key, value in text_batch.items()})
    image_loader = DataLoader(ImageDataset(train, image_transform()), batch_size=4, shuffle=False, num_workers=0)
    image_model = create_resnet().to(device)
    image_batch = next(iter(image_loader))
    with torch.no_grad(), torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
        image_logits = image_model(image_batch["image"].to(device))
    if text_out.logits.shape != (8, 2) or image_logits.shape != (4, 2):
        raise ValueError("Unexpected smoke-test output shape")
    if not np.array_equal(text_batch["labels"].numpy(), train.iloc[text_indices.numpy()]["label"].to_numpy()):
        raise ValueError("Text labels are not aligned")
    if not np.array_equal(image_batch["label"].numpy(), train.iloc[image_batch["sample_index"].numpy()]["label"].to_numpy()):
        raise ValueError("Image labels are not aligned")
    result = {"passed": True, "device": str(device), "gpu": torch.cuda.get_device_name(0) if device.type == "cuda" else None, "text_batch_shape": list(text_out.logits.shape), "image_batch_shape": list(image_logits.shape), "labels_aligned": True, "output_root": str(root)}
    dump_json(paths(root)["logs"] / "smoke_test.json", result)
    print(json.dumps(result, indent=2))


def train_roberta(root: Path, epochs: int, batch_size: int) -> None:
    p = paths(root)
    if (p["roberta_checkpoint"] / "model.safetensors").exists() or (p["roberta_checkpoint"] / "pytorch_model.bin").exists():
        raise FileExistsError("RoBERTa checkpoint already exists; refusing to overwrite it")
    set_seed()
    df = load_manifest(root)
    train, validation = split_df(df, "train"), split_df(df, "validation")
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    tokenizer = AutoTokenizer.from_pretrained(MODEL_NAME)
    train_loader = DataLoader(TextDataset(train, tokenizer), batch_size=batch_size, shuffle=True, num_workers=0, pin_memory=device.type == "cuda", generator=torch.Generator().manual_seed(SEED))
    validation_loader = DataLoader(TextDataset(validation, tokenizer), batch_size=batch_size, shuffle=False, num_workers=0, pin_memory=device.type == "cuda")
    model = AutoModelForSequenceClassification.from_pretrained(MODEL_NAME, num_labels=2).to(device)
    optimizer = AdamW(model.parameters(), lr=2e-5, weight_decay=0.01)
    total_steps = len(train_loader) * epochs
    scheduler = get_linear_schedule_with_warmup(optimizer, num_warmup_steps=int(total_steps * 0.10), num_training_steps=total_steps)
    scaler = torch.amp.GradScaler("cuda", enabled=device.type == "cuda")
    history, best = [], -1.0
    for epoch in range(1, epochs + 1):
        model.train()
        total_loss = 0.0
        for step, batch in enumerate(train_loader, 1):
            batch.pop("sample_index")
            batch = {key: value.to(device, non_blocking=True) for key, value in batch.items()}
            optimizer.zero_grad(set_to_none=True)
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                output = model(**batch)
                loss = output.loss
            scaler.scale(loss).backward()
            scaler.unscale_(optimizer)
            torch.nn.utils.clip_grad_norm_(model.parameters(), 1.0)
            scaler.step(optimizer)
            scaler.update()
            scheduler.step()
            total_loss += float(loss.item())
            if step % 100 == 0:
                print(f"RoBERTa epoch {epoch} step {step}/{len(train_loader)} loss={total_loss/step:.4f}", flush=True)
        val_metrics, indices, labels, preds, probs = text_evaluate(model, validation_loader, device)
        record = {"epoch": epoch, "train_loss": total_loss / len(train_loader), **{f"validation_{k}": v for k, v in val_metrics.items() if k != "confusion_matrix"}}
        history.append(record)
        print(json.dumps(record, allow_nan=False), flush=True)
        if val_metrics["macro_f1"] > best:
            best = val_metrics["macro_f1"]
            model.save_pretrained(p["roberta_checkpoint"])
            tokenizer.save_pretrained(p["roberta_checkpoint"])
            prediction_frame(validation, indices, labels, preds, probs, "roberta").to_csv(p["predictions"] / "roberta_validation.csv", index=False)
            dump_json(p["metrics"] / "roberta_best_validation.json", {"best_epoch": epoch, "metrics": val_metrics, "checkpoint": str(p["roberta_checkpoint"])})
    pd.DataFrame(history).to_csv(p["metrics"] / "roberta_training_history.csv", index=False)
    print(f"Best validation macro F1: {best:.6f}")


def train_resnet(root: Path, epochs: int, batch_size: int, num_workers: int) -> None:
    p = paths(root)
    checkpoint_path = p["resnet_checkpoint"] / "best_model.pt"
    if checkpoint_path.exists():
        raise FileExistsError("ResNet checkpoint already exists; refusing to overwrite it")
    set_seed()
    df = load_manifest(root)
    train, validation = split_df(df, "train"), split_df(df, "validation")
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    loader_args = {"num_workers": num_workers, "pin_memory": device.type == "cuda", "worker_init_fn": worker_seed}
    if num_workers > 0:
        loader_args["persistent_workers"] = True
    train_loader = DataLoader(ImageDataset(train, image_transform()), batch_size=batch_size, shuffle=True, generator=torch.Generator().manual_seed(SEED), **loader_args)
    validation_loader = DataLoader(ImageDataset(validation, image_transform()), batch_size=batch_size, shuffle=False, **loader_args)
    model = create_resnet().to(device)
    criterion = nn.CrossEntropyLoss()
    optimizer = AdamW(model.parameters(), lr=1e-4, weight_decay=0.01)
    scaler = torch.amp.GradScaler("cuda", enabled=device.type == "cuda")
    history, best = [], -1.0
    for epoch in range(1, epochs + 1):
        model.train()
        total_loss = 0.0
        for step, batch in enumerate(train_loader, 1):
            images = batch["image"].to(device, non_blocking=True)
            labels = batch["label"].to(device, non_blocking=True)
            optimizer.zero_grad(set_to_none=True)
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                logits = model(images)
                loss = criterion(logits, labels)
            scaler.scale(loss).backward()
            scaler.unscale_(optimizer)
            torch.nn.utils.clip_grad_norm_(model.parameters(), 1.0)
            scaler.step(optimizer)
            scaler.update()
            total_loss += float(loss.item())
            if step % 50 == 0:
                print(f"ResNet epoch {epoch} step {step}/{len(train_loader)} loss={total_loss/step:.4f}", flush=True)
        val_metrics, indices, labels, preds, probs = image_evaluate(model, validation_loader, device)
        record = {"epoch": epoch, "train_loss": total_loss / len(train_loader), **{f"validation_{k}": v for k, v in val_metrics.items() if k != "confusion_matrix"}}
        history.append(record)
        print(json.dumps(record, allow_nan=False), flush=True)
        if val_metrics["macro_f1"] > best:
            best = val_metrics["macro_f1"]
            torch.save({"model_state_dict": model.state_dict(), "model": "resnet50", "weights": "IMAGENET1K_V2", "num_classes": 2, "best_epoch": epoch, "validation_macro_f1": best}, checkpoint_path)
            prediction_frame(validation, indices, labels, preds, probs, "resnet").to_csv(p["predictions"] / "resnet_validation.csv", index=False)
            dump_json(p["metrics"] / "resnet_best_validation.json", {"best_epoch": epoch, "metrics": val_metrics, "checkpoint": str(checkpoint_path)})
    pd.DataFrame(history).to_csv(p["metrics"] / "resnet_training_history.csv", index=False)
    print(f"Best validation macro F1: {best:.6f}")


def stage_lock(root: Path) -> None:
    p = paths(root)
    if p["lock"].exists():
        raise FileExistsError("Validation lock already exists; refusing to replace it")
    text = pd.read_csv(p["predictions"] / "roberta_validation.csv")
    image = pd.read_csv(p["predictions"] / "resnet_validation.csv")
    merged = text.merge(image, on=["sample_id", "true_label"], validate="one_to_one")
    expected = len(split_df(load_manifest(root), "validation"))
    if len(merged) != expected:
        raise ValueError(f"Paired validation count {len(merged)} does not equal {expected}")
    merged.to_csv(p["predictions"] / "validation_predictions.csv", index=False)
    rows = []
    y = merged["true_label"].to_numpy(dtype=int)
    for alpha in np.arange(0, 1.0001, 0.05):
        probability = alpha * merged["roberta_probability_class1"].to_numpy() + (1 - alpha) * merged["resnet_probability_class1"].to_numpy()
        pred = (probability >= THRESHOLD).astype(int)
        score = metrics_for(y, pred, probability)
        rows.append({"alpha_text": round(float(alpha), 2), "alpha_image": round(float(1-alpha), 2), **{k: v for k, v in score.items() if k not in {"confusion_matrix", "recall_class_0", "recall_class_1"}}})
    search = pd.DataFrame(rows)
    search.to_csv(p["metrics"] / "validation_alpha_search.csv", index=False)
    maximum = search["macro_f1"].max()
    tied = search[np.isclose(search["macro_f1"], maximum)].copy()
    tied["distance_from_half"] = (tied["alpha_text"] - 0.5).abs()
    selected = tied.sort_values(["distance_from_half", "alpha_text"], ascending=[True, True]).iloc[0]

    # Optional fair text control: tune threshold and Platt calibration on validation only.
    threshold_rows = []
    for threshold in np.arange(0.05, 0.951, 0.01):
        pred = (merged["roberta_probability_class1"].to_numpy() >= threshold).astype(int)
        threshold_rows.append({"threshold": round(float(threshold), 2), "macro_f1": f1_score(y, pred, average="macro", zero_division=0)})
    threshold_search = pd.DataFrame(threshold_rows)
    threshold_search.to_csv(p["metrics"] / "roberta_validation_threshold_search.csv", index=False)
    threshold_best = threshold_search.sort_values(["macro_f1", "threshold"], ascending=[False, True]).iloc[0]
    calibrator = LogisticRegression(random_state=SEED).fit(merged[["roberta_probability_class1"]], y)
    dump_json(p["metrics"] / "fair_text_validation_control.json", {"selected_threshold": float(threshold_best["threshold"]), "validation_macro_f1": float(threshold_best["macro_f1"]), "platt_coefficient": float(calibrator.coef_[0, 0]), "platt_intercept": float(calibrator.intercept_[0])})

    lock = {"locked_utc": datetime.now(timezone.utc).isoformat(), "selection_partition": "validation", "paired_validation_samples": int(len(merged)), "selection_metric": "macro_f1", "selected_alpha_text": float(selected["alpha_text"]), "selected_alpha_image": float(selected["alpha_image"]), "validation_macro_f1": float(selected["macro_f1"]), "classification_threshold": THRESHOLD, "tied_alpha_values": tied["alpha_text"].astype(float).tolist(), "tie_break": "closest to 0.50, then lower alpha", "roberta_checkpoint": str(p["roberta_checkpoint"]), "resnet_checkpoint": str(p["resnet_checkpoint"] / "best_model.pt")}
    dump_json(p["lock"], lock)
    config = json.loads(p["config"].read_text(encoding="utf-8"))
    config["fusion"]["selected_alpha"] = lock["selected_alpha_text"]
    config["fusion"]["locked_utc"] = lock["locked_utc"]
    dump_json(p["config"], config)
    print(json.dumps(lock, indent=2))


# END REGISTERED SOURCE BLOCK


In [88]:
%%project_source v2/experiments/source_disjoint/run_source_disjoint.py 3
def ece(labels, probabilities, n_bins=N_BINS):
    labels = np.asarray(labels, dtype=int)
    probabilities = np.asarray(probabilities, dtype=float)
    predictions = (probabilities >= 0.5).astype(int)
    confidence = np.maximum(probabilities, 1 - probabilities)
    correctness = (predictions == labels).astype(float)
    edges = np.linspace(0.5, 1.0, n_bins + 1)
    value, rows = 0.0, []
    for index, (lower, upper) in enumerate(zip(edges[:-1], edges[1:])):
        mask = (confidence >= lower) & (confidence <= upper if index == n_bins - 1 else confidence < upper)
        count = int(mask.sum())
        mean_confidence = float(confidence[mask].mean()) if count else None
        accuracy = float(correctness[mask].mean()) if count else None
        gap = abs(accuracy - mean_confidence) if count else None
        if count:
            value += count / len(labels) * gap
        rows.append({"bin_lower": float(lower), "bin_upper": float(upper), "count": count, "mean_confidence": mean_confidence, "accuracy": accuracy, "gap": gap})
    return float(value), rows


def calibration_for(name, labels, probabilities):
    clipped = np.clip(np.asarray(probabilities, dtype=float), 1e-7, 1 - 1e-7)
    ece_value, bins = ece(labels, clipped)
    return {"model": name, "brier": float(brier_score_loss(labels, clipped)), "log_loss": float(log_loss(labels, clipped)), "ece": ece_value}, bins


def bootstrap(root: Path, y, models: dict[str, tuple[np.ndarray, np.ndarray]]) -> pd.DataFrame:
    rng = np.random.default_rng(SEED)
    text_pred, text_prob = models["roberta"]
    fusion_pred, fusion_prob = models["late_fusion"]
    observed_text = metrics_for(y, text_pred, text_prob)
    observed_fusion = metrics_for(y, fusion_pred, fusion_prob)
    names = ["accuracy", "f1", "macro_f1", "roc_auc", "pr_auc"]
    values = {name: [] for name in names}
    for _ in range(N_BOOTSTRAPS):
        idx = rng.integers(0, len(y), size=len(y))
        ys = y[idx]
        basic_text = metrics_for(ys, text_pred[idx], text_prob[idx])
        basic_fusion = metrics_for(ys, fusion_pred[idx], fusion_prob[idx])
        for name in names:
            if basic_text[name] is not None and basic_fusion[name] is not None:
                values[name].append(basic_fusion[name] - basic_text[name])
    pd.DataFrame({name: pd.Series(series) for name, series in values.items()}).to_csv(paths(root)["bootstrap"] / "paired_differences.csv", index=False)
    rows = []
    for name in names:
        series = np.asarray(values[name])
        rows.append({"metric": name, "difference": observed_fusion[name] - observed_text[name], "ci_lower": float(np.percentile(series, 2.5)), "ci_upper": float(np.percentile(series, 97.5)), "valid_iterations": int(len(series)), "requested_iterations": N_BOOTSTRAPS})
    result = pd.DataFrame(rows)
    result.to_csv(paths(root)["metrics"] / "statistical_comparison.csv", index=False)
    return result


def reliability_plot(root: Path, bins_by_model: dict[str, list[dict]]) -> None:
    fig, ax = plt.subplots(figsize=(7, 6))
    ax.plot([0.5, 1.0], [0.5, 1.0], color="black", linestyle=":", label="Perfect calibration")
    for name, rows in bins_by_model.items():
        frame = pd.DataFrame(rows).dropna(subset=["mean_confidence", "accuracy"])
        ax.plot(frame["mean_confidence"], frame["accuracy"], marker="o", label=name)
    ax.set(xlabel="Mean confidence", ylabel="Observed accuracy", xlim=(0.5, 1.0), ylim=(0.5, 1.0), title="Source-disjoint test reliability")
    ax.legend()
    fig.tight_layout()
    fig.savefig(paths(root)["figures"] / "reliability_diagram.png", dpi=180)
    plt.close(fig)


def markdown_table(frame: pd.DataFrame, decimals: int = 4) -> str:
    """Render a small DataFrame without the optional tabulate dependency."""
    display = frame.copy()
    for column in display.select_dtypes(include=["float", "floating"]).columns:
        display[column] = display[column].map(lambda value: "" if pd.isna(value) else f"{value:.{decimals}f}")
    headers = [str(column) for column in display.columns]
    lines = ["| " + " | ".join(headers) + " |", "| " + " | ".join(["---"] * len(headers)) + " |"]
    for row in display.itertuples(index=False, name=None):
        lines.append("| " + " | ".join(str(value).replace("|", "\\|") for value in row) + " |")
    return "\n".join(lines)


def stage_test(root: Path, text_batch: int, image_batch: int, num_workers: int) -> None:
    p = paths(root)
    final_predictions_path = p["predictions"] / "test_predictions.csv"
    if final_predictions_path.exists():
        raise FileExistsError("Test predictions already exist; refusing to evaluate the locked test twice")
    lock = json.loads(p["lock"].read_text(encoding="utf-8"))
    alpha = float(lock["selected_alpha_text"])
    set_seed()
    test = split_df(load_manifest(root), "test")
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")

    tokenizer = AutoTokenizer.from_pretrained(p["roberta_checkpoint"])
    text_loader = DataLoader(TextDataset(test, tokenizer), batch_size=text_batch, shuffle=False, num_workers=0, pin_memory=device.type == "cuda")
    text_model = AutoModelForSequenceClassification.from_pretrained(p["roberta_checkpoint"]).to(device)
    _, ti, ty, tp, tprob = text_evaluate(text_model, text_loader, device)
    text_frame = prediction_frame(test, ti, ty, tp, tprob, "roberta")
    del text_model
    if device.type == "cuda":
        torch.cuda.empty_cache()

    loader_args = {"num_workers": num_workers, "pin_memory": device.type == "cuda", "worker_init_fn": worker_seed}
    if num_workers > 0:
        loader_args["persistent_workers"] = True
    image_loader = DataLoader(ImageDataset(test, image_transform()), batch_size=image_batch, shuffle=False, **loader_args)
    image_model = create_resnet().to(device)
    checkpoint = torch.load(p["resnet_checkpoint"] / "best_model.pt", map_location=device, weights_only=True)
    image_model.load_state_dict(checkpoint["model_state_dict"])
    _, ii, iy, ip, iprob = image_evaluate(image_model, image_loader, device)
    image_frame = prediction_frame(test, ii, iy, ip, iprob, "resnet")

    predictions = text_frame.merge(image_frame, on=["sample_id", "true_label"], validate="one_to_one")
    diagnostics = test[["id", "subreddit"]].rename(columns={"id": "sample_id"})
    predictions = predictions.merge(diagnostics, on="sample_id", validate="one_to_one")
    predictions["fusion_probability_class1"] = alpha * predictions["roberta_probability_class1"] + (1 - alpha) * predictions["resnet_probability_class1"]
    predictions["fusion_prediction"] = (predictions["fusion_probability_class1"] >= THRESHOLD).astype(int)
    predictions.to_csv(final_predictions_path, index=False)

    y = predictions["true_label"].to_numpy(dtype=int)
    model_arrays = {
        "roberta": (predictions["roberta_prediction"].to_numpy(dtype=int), predictions["roberta_probability_class1"].to_numpy()),
        "resnet50": (predictions["resnet_prediction"].to_numpy(dtype=int), predictions["resnet_probability_class1"].to_numpy()),
        "late_fusion": (predictions["fusion_prediction"].to_numpy(dtype=int), predictions["fusion_probability_class1"].to_numpy()),
    }
    metric_rows, full_metrics = [], {}
    calibration_rows, bins_by_model = [], {}
    for name, (pred, prob) in model_arrays.items():
        values = metrics_for(y, pred, prob)
        full_metrics[name] = values
        cal, bins = calibration_for(name, y, prob)
        calibration_rows.append(cal)
        bins_by_model[name] = bins
        pd.DataFrame(bins).to_csv(p["calibration"] / f"{name}_bins.csv", index=False)
        metric_rows.append({"model": name, **{key: value for key, value in values.items() if key != "confusion_matrix"}, **{key: value for key, value in cal.items() if key != "model"}})
    metric_summary = pd.DataFrame(metric_rows)
    metric_summary.to_csv(p["metrics"] / "summary.csv", index=False)
    dump_json(p["metrics"] / "summary.json", {"test_samples": len(predictions), "selected_alpha_text": alpha, "models": full_metrics})
    calibration_frame = pd.DataFrame(calibration_rows)
    calibration_frame.to_csv(p["calibration"] / "calibration_metrics.csv", index=False)
    dump_json(p["calibration"] / "calibration_metrics.json", {"n_bins": N_BINS, "convention": "confidence bins from 0.5 to 1.0", "models": calibration_rows})
    reliability_plot(root, bins_by_model)

    cr = model_arrays["roberta"][0] == y
    ci = model_arrays["resnet50"][0] == y
    cf = model_arrays["late_fusion"][0] == y
    b = int(np.sum(cr & ~cf))
    c = int(np.sum(~cr & cf))
    mcnemar_p = float(binomtest(min(b, c), n=b + c, p=0.5, alternative="two-sided").pvalue) if b + c else 1.0
    mcnemar = {"both_correct": int(np.sum(cr & cf)), "both_wrong": int(np.sum(~cr & ~cf)), "roberta_correct_fusion_wrong": b, "fusion_correct_roberta_wrong": c, "discordant": b + c, "exact_p_value": mcnemar_p}
    dump_json(p["metrics"] / "mcnemar.json", mcnemar)
    stats = bootstrap(root, y, model_arrays)
    complementarity = {
        "roberta_vs_fusion": mcnemar,
        "roberta_vs_resnet_disagreements": int(np.sum(model_arrays["roberta"][0] != model_arrays["resnet50"][0])),
        "roberta_only_correct": int(np.sum(cr & ~ci)),
        "resnet_only_correct": int(np.sum(~cr & ci)),
        "image_correct_text_wrong_recovered_by_fusion": int(np.sum(~cr & ci & cf)),
        "text_correct_image_wrong_preserved_by_fusion": int(np.sum(cr & ~ci & cf)),
    }
    dump_json(p["metrics"] / "error_complementarity.json", complementarity)

    # Apply the validation-selected fair text threshold and Platt model once to test.
    fair = json.loads((p["metrics"] / "fair_text_validation_control.json").read_text(encoding="utf-8"))
    tuned_pred = (model_arrays["roberta"][1] >= fair["selected_threshold"]).astype(int)
    z = fair["platt_intercept"] + fair["platt_coefficient"] * model_arrays["roberta"][1]
    platt_prob = 1 / (1 + np.exp(-z))
    pd.DataFrame([
        {"control": "validation_tuned_threshold", "threshold": fair["selected_threshold"], **{k: v for k, v in metrics_for(y, tuned_pred, model_arrays["roberta"][1]).items() if k != "confusion_matrix"}},
        {"control": "validation_platt_calibration", "threshold": 0.5, **{k: v for k, v in metrics_for(y, (platt_prob >= 0.5).astype(int), platt_prob).items() if k != "confusion_matrix"}},
    ]).to_csv(p["metrics"] / "fair_text_test_control.csv", index=False)

    original = {"roberta": {"accuracy": 0.8046, "macro_f1": 0.8000, "roc_auc": 0.8846, "pr_auc": 0.9027}, "resnet50": {"accuracy": 0.7382, "macro_f1": 0.7275, "roc_auc": 0.7976, "pr_auc": 0.8053}, "late_fusion": {"accuracy": 0.8242, "macro_f1": 0.8188, "roc_auc": 0.8993, "pr_auc": 0.9097}}
    penalty_rows = []
    for name in original:
        for metric, old in original[name].items():
            penalty_rows.append({"model": name, "metric": metric, "ordinary_locked_holdout": old, "source_disjoint": full_metrics[name][metric], "change_source_disjoint_minus_ordinary": full_metrics[name][metric] - old})
    pd.DataFrame(penalty_rows).to_csv(p["metrics"] / "generalisation_penalty.csv", index=False)

    counts = pd.read_csv(p["manifests"] / "split_counts.csv")
    macro_row = stats[stats["metric"].eq("macro_f1")].iloc[0]
    best_text = json.loads((p["metrics"] / "roberta_best_validation.json").read_text(encoding="utf-8"))
    best_image = json.loads((p["metrics"] / "resnet_best_validation.json").read_text(encoding="utf-8"))
    lines = [
        "# Source-disjoint evaluation results", "",
        "## Dataset and split verification", "",
        "The manifest assigns every subreddit to one partition. No subreddit appears in more than one split. Both labels occur in every split. All image files opened correctly and the known regional-unavailable placeholder was absent.", "",
        markdown_table(counts), "",
        "The source-disjoint manifest was created from the existing cleaned multimodal pool. The manifest count is therefore also the final usable count, with no further removals in this run.", "",
        "## Locked validation choices", "",
        f"RoBERTa checkpoint: `{best_text['checkpoint']}` (epoch {best_text['best_epoch']}).", "",
        f"ResNet-50 checkpoint: `{best_image['checkpoint']}` (epoch {best_image['best_epoch']}).", "",
        f"Validation selected alpha = {alpha:.2f} for RoBERTa and {1-alpha:.2f} for ResNet-50. The classification threshold remained 0.50.", "",
        "The complete search is in `metrics/validation_alpha_search.csv`.", "",
        "## Source-disjoint test performance", "", markdown_table(metric_summary), "",
        "## Calibration", "", markdown_table(calibration_frame), "",
        "Lower Brier score, log loss and ECE indicate better calibration.", "",
        "## Paired statistical comparison", "",
        f"Late fusion and RoBERTa were compared on {len(y):,} paired test cases. Both were correct on {mcnemar['both_correct']:,}; both were wrong on {mcnemar['both_wrong']:,}. RoBERTa alone was correct on {b:,} and fusion alone on {c:,}. The exact McNemar p-value was {mcnemar_p:.6g}.", "",
        markdown_table(stats), "",
        "## Error complementarity", "",
        f"RoBERTa and ResNet-50 disagreed on {complementarity['roberta_vs_resnet_disagreements']:,} cases. RoBERTa alone was correct on {complementarity['roberta_only_correct']:,}; ResNet-50 alone was correct on {complementarity['resnet_only_correct']:,}. Late fusion recovered {complementarity['image_correct_text_wrong_recovered_by_fusion']:,} image-correct/text-wrong cases and preserved {complementarity['text_correct_image_wrong_preserved_by_fusion']:,} text-correct/image-wrong cases.", "",
        "## Interpretation", "",
        f"Removing subreddit overlap changed RoBERTa macro F1 by {full_metrics['roberta']['macro_f1']-0.8000:+.4f}, ResNet-50 by {full_metrics['resnet50']['macro_f1']-0.7275:+.4f}, and late fusion by {full_metrics['late_fusion']['macro_f1']-0.8188:+.4f} compared with the ordinary locked holdout. Late fusion changed macro F1 over RoBERTa by {full_metrics['late_fusion']['macro_f1']-full_metrics['roberta']['macro_f1']:+.4f}. Its paired 95% bootstrap interval was [{macro_row['ci_lower']:+.4f}, {macro_row['ci_upper']:+.4f}]. Validation selected zero text weight, so the locked late-fusion result is identical to ResNet-50 and does not show a benefit from combining modalities. These figures measure transfer to unseen subreddit groups rather than performance on the earlier mixed-source holdout.", "",
    ]
    (p["reports"] / "source_disjoint_results.md").write_text("\n".join(lines), encoding="utf-8")
    config = json.loads(p["config"].read_text(encoding="utf-8"))
    config["test_evaluated_utc"] = datetime.now(timezone.utc).isoformat()
    config["test_predictions"] = str(final_predictions_path)
    dump_json(p["config"], config)
    print(metric_summary.to_string(index=False))
    print(json.dumps(mcnemar, indent=2))


# END REGISTERED SOURCE BLOCK


In [89]:
%%project_source v2/experiments/source_disjoint/run_source_disjoint.py 4
def main() -> None:
    parser = argparse.ArgumentParser()
    parser.add_argument("stage", choices=["audit", "smoke", "train-roberta", "train-resnet", "lock", "test"])
    parser.add_argument("--experiment-root", type=Path, default=DEFAULT_EXPERIMENT_ROOT)
    parser.add_argument("--epochs", type=int, default=3)
    parser.add_argument("--batch-size", type=int)
    parser.add_argument("--num-workers", type=int, default=2)
    args = parser.parse_args()
    root = args.experiment_root.resolve()
    if args.stage == "audit": stage_audit(root)
    elif args.stage == "smoke": stage_smoke(root)
    elif args.stage == "train-roberta": train_roberta(root, args.epochs, args.batch_size or 16)
    elif args.stage == "train-resnet": train_resnet(root, args.epochs, args.batch_size or 32, args.num_workers)
    elif args.stage == "lock": stage_lock(root)
    elif args.stage == "test": stage_test(root, args.batch_size or 16, 32, args.num_workers)


if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


<a id="support"></a>
## 10. Verification, configuration and historical sources

### 10.1 Verify saved results

Verify archived evidence fingerprints and recompute headline metrics from saved predictions without running model inference.

**Source:** `tools/verify_saved_results.py`  
**Imported modules:** `csv`, `hashlib`, `json`, `math`, `pathlib`  
**Top-level components:** `require`, `load_csv`, `verify_models`, `main`

The following cells contain the complete source; Run All registers it for inspection/export.

In [90]:
%%project_source tools/verify_saved_results.py 0
"""Read-only verification of the packaged dissertation evidence (stdlib only)."""
from pathlib import Path
import csv
import hashlib
import json
import math

ROOT = Path(__file__).resolve().parents[1]


def require(condition, message):
    if not condition:
        raise AssertionError(message)


def load_csv(path):
    with path.open(encoding="utf-8-sig", newline="") as handle:
        return list(csv.DictReader(handle))


def verify_models(rows, label, specs, scores, macro_key):
    for model, prediction, probability in specs:
        cm = [[0, 0], [0, 0]]
        for row in rows:
            y, pred, prob = int(row[label]), int(row[prediction]), float(row[probability])
            require(y in (0, 1) and pred in (0, 1), "Invalid binary label")
            require(math.isfinite(prob) and 0 <= prob <= 1, "Invalid probability")
            require(pred == int(prob >= 0.5), f"{model}: prediction/threshold mismatch")
            cm[y][pred] += 1
        accuracy = (cm[0][0] + cm[1][1]) / len(rows)
        macro = sum(2 * cm[k][k] / (2 * cm[k][k] + cm[0][1] + cm[1][0]) for k in (0, 1)) / 2
        require(cm == scores[model]["confusion_matrix"], f"{model}: confusion matrix mismatch")
        require(abs(accuracy - scores[model]["accuracy"]) < 1e-10, f"{model}: accuracy mismatch")
        require(abs(macro - scores[model][macro_key]) < 1e-10, f"{model}: macro F1 mismatch")
        print(f"  {model:12s} n={len(rows):4d} accuracy={accuracy:.4f} macro_F1={macro:.4f}")


def main():
    manifest = load_csv(ROOT / "evidence_manifest.csv")
    for row in manifest:
        path = ROOT / row["path"]
        require(path.is_file(), f"Missing evidence: {row['path']}")
        require(path.stat().st_size == int(row["bytes"]), f"Size changed: {row['path']}")
        require(hashlib.sha256(path.read_bytes()).hexdigest() == row["sha256"], f"Fingerprint changed: {row['path']}")
    print(f"Verified {len(manifest)} evidence fingerprints.")

    ordinary = ROOT / "multimodal-fake-news-detection/results/metrics/final_evaluation"
    rows = load_csv(ordinary / "final_predictions.csv")
    saved = json.loads((ordinary / "final_results.json").read_text())
    ids = [r["id"] for r in rows]
    require(len(ids) == len(set(ids)) == saved["holdout"]["samples"] == 5000, "Ordinary ID/size mismatch")
    require(hashlib.sha256("\n".join(ids).encode()).hexdigest() == saved["holdout"]["ordered_id_sha256"], "Ordinary ordered-ID freeze mismatch")
    alpha = saved["locked_specification"]["alpha_text"]
    require(alpha == 0.45, "Unexpected ordinary fusion weight")
    for r in rows:
        expected = alpha * float(r["probability_roberta"]) + (1-alpha) * float(r["probability_resnet"])
        require(abs(expected-float(r["probability_fusion"])) < 1e-10, "Ordinary fusion arithmetic mismatch")
    print("Ordinary locked holdout:")
    verify_models(rows, "label", [(m, f"prediction_{col}", f"probability_{col}") for m,col in [("roberta","roberta"),("resnet","resnet"),("late_fusion","fusion")]], saved["metrics"], "f1_macro")

    source = ROOT / "v2/experiments/source_disjoint"
    rows = load_csv(source / "predictions/test_predictions.csv")
    saved = json.loads((source / "metrics/summary.json").read_text())
    require(len(rows) == len({r["sample_id"] for r in rows}) == saved["test_samples"] == 2739, "Source ID/size mismatch")
    require(saved["selected_alpha_text"] == 0, "Unexpected source-disjoint weight")
    for r in rows:
        require(abs(float(r["fusion_probability_class1"])-float(r["resnet_probability_class1"])) < 1e-10, "Source fusion arithmetic mismatch")
    print("Source-disjoint test:")
    verify_models(rows, "true_label", [(m, f"{col}_prediction", f"{col}_probability_class1") for m,col in [("roberta","roberta"),("resnet50","resnet"),("late_fusion","fusion")]], saved["models"], "macro_f1")
    print("PASS: packaged results agree with saved predictions. No experiments were rerun.")


if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


### 10.2 Test environment

Project support implementation.

**Source:** `multimodal-fake-news-detection/tests/test_environment.py`  
**Imported modules:** `torch`  
**Top-level components:** `test_pytorch_available`, `test_tensor_creation`

The following cells contain the complete source; Run All registers it for inspection/export.

In [91]:
%%project_source multimodal-fake-news-detection/tests/test_environment.py 0
import torch


def test_pytorch_available():
    assert torch.__version__ is not None


def test_tensor_creation():
    tensor = torch.tensor([1.0, 2.0, 3.0])
    assert tensor.shape == (3,)
# END REGISTERED SOURCE BLOCK


### Package module: `multimodal-fake-news-detection/src/fake_news/__init__.py`

Preserved even where it is an empty package initialiser.

In [92]:
%%project_source multimodal-fake-news-detection/src/fake_news/__init__.py 0

# END REGISTERED SOURCE BLOCK


### Package module: `multimodal-fake-news-detection/src/fake_news/data/__init__.py`

Preserved even where it is an empty package initialiser.

In [93]:
%%project_source multimodal-fake-news-detection/src/fake_news/data/__init__.py 0

# END REGISTERED SOURCE BLOCK


### Package module: `multimodal-fake-news-detection/src/fake_news/evaluation/__init__.py`

Preserved even where it is an empty package initialiser.

In [94]:
%%project_source multimodal-fake-news-detection/src/fake_news/evaluation/__init__.py 0

# END REGISTERED SOURCE BLOCK


### Package module: `multimodal-fake-news-detection/src/fake_news/explainability/__init__.py`

Preserved even where it is an empty package initialiser.

In [95]:
%%project_source multimodal-fake-news-detection/src/fake_news/explainability/__init__.py 0

# END REGISTERED SOURCE BLOCK


### Package module: `multimodal-fake-news-detection/src/fake_news/models/__init__.py`

Preserved even where it is an empty package initialiser.

In [96]:
%%project_source multimodal-fake-news-detection/src/fake_news/models/__init__.py 0

# END REGISTERED SOURCE BLOCK


### Package module: `multimodal-fake-news-detection/src/fake_news/training/__init__.py`

Preserved even where it is an empty package initialiser.

In [97]:
%%project_source multimodal-fake-news-detection/src/fake_news/training/__init__.py 0

# END REGISTERED SOURCE BLOCK


### Historical local variants

These are provenance copies, not extra experiments. The local source-disjoint runner and report builder contain hard-coded F: paths; the runner helper below refuses to execute anything under `historical/`. Use the canonical runner for reproduction. The earlier methodology setup is also retained. Other local Python scripts were compared with the submission copy and were identical.

#### Earlier local file: `v2/experiments/source_disjoint/run_source_disjoint.py`

In [98]:
%%project_source historical/v2/experiments/source_disjoint/run_source_disjoint.py 0
"""Isolated source-disjoint retraining and evaluation for the Fakeddit study.

The command is deliberately split into stages so the test partition is not used
until both validation checkpoints and the late-fusion coefficient are locked.
"""

from __future__ import annotations

import argparse
import hashlib
import json
import os
import platform
import random
import shutil
import sys
from datetime import datetime, timezone
from pathlib import Path

import matplotlib.pyplot as plt
import numpy as np
import pandas as pd
import scipy
import sklearn
import torch
import torch.nn as nn
import torchvision
import transformers
from PIL import Image
from scipy.stats import binomtest
from sklearn.linear_model import LogisticRegression
from sklearn.metrics import (
    accuracy_score,
    average_precision_score,
    brier_score_loss,
    confusion_matrix,
    f1_score,
    log_loss,
    precision_score,
    recall_score,
    roc_auc_score,
)
from torch.optim import AdamW
from torch.utils.data import DataLoader, Dataset
from torchvision import transforms
from torchvision.models import ResNet50_Weights, resnet50
from transformers import (
    AutoModelForSequenceClassification,
    AutoTokenizer,
    get_linear_schedule_with_warmup,
)


SEED = 42
MODEL_NAME = "roberta-base"
MAX_LENGTH = 64
THRESHOLD = 0.50
N_BINS = 10
N_BOOTSTRAPS = 5000
PLACEHOLDER_SHA256 = "faa24ec881e6040655c187a681d6dc496eb8aa41e1bd0652a180b3a40b457187"
PROJECT_ROOT = Path(r"F:\data sci\project\multimodal-fake-news-detection")
SOURCE_MANIFEST = Path(r"F:\data sci\project\v2\manifests\source_disjoint.parquet")
DEFAULT_EXPERIMENT_ROOT = Path(r"F:\data sci\project\v2\experiments\source_disjoint")


def paths(root: Path) -> dict[str, Path]:
    return {
        "root": root,
        "manifests": root / "manifests",
        "checkpoints": root / "checkpoints",
        "roberta_checkpoint": root / "checkpoints" / "roberta",
        "resnet_checkpoint": root / "checkpoints" / "resnet50",
        "predictions": root / "predictions",
        "metrics": root / "metrics",
        "logs": root / "logs",
        "figures": root / "figures",
        "bootstrap": root / "bootstrap",
        "calibration": root / "calibration",
        "reports": root / "reports",
        "manifest": root / "manifests" / "source_disjoint.parquet",
        "config": root / "experiment_config.json",
        "audit": root / "manifests" / "manifest_audit.json",
        "lock": root / "metrics" / "validation_lock.json",
    }


def make_dirs(root: Path) -> None:
    for key, value in paths(root).items():
        if key not in {"manifest", "config", "audit", "lock"}:
            value.mkdir(parents=True, exist_ok=True)


def dump_json(path: Path, value: dict) -> None:
    path.parent.mkdir(parents=True, exist_ok=True)
    path.write_text(json.dumps(value, indent=2, allow_nan=False), encoding="utf-8")


def set_seed(seed: int = SEED) -> None:
    os.environ["PYTHONHASHSEED"] = str(seed)
    random.seed(seed)
    np.random.seed(seed)
    torch.manual_seed(seed)
    if torch.cuda.is_available():
        torch.cuda.manual_seed_all(seed)
    torch.backends.cudnn.deterministic = True
    torch.backends.cudnn.benchmark = False


def resolve_image_path(value: str) -> Path:
    path = Path(str(value))
    return path if path.is_absolute() else PROJECT_ROOT / path


def load_manifest(root: Path) -> pd.DataFrame:
    path = paths(root)["manifest"]
    if not path.exists():
        raise FileNotFoundError(f"Run the audit stage first: {path}")
    df = pd.read_parquet(path)
    required = {"id", "label", "text", "image_path", "subreddit", "v2_split"}
    missing = required.difference(df.columns)
    if missing:
        raise ValueError(f"Manifest lacks columns: {sorted(missing)}")
    df = df.copy()
    df["id"] = df["id"].astype(str)
    df["label"] = df["label"].astype(int)
    df["resolved_image_path"] = df["image_path"].map(lambda x: str(resolve_image_path(x)))
    return df


def split_df(df: pd.DataFrame, split: str) -> pd.DataFrame:
    result = df.loc[df["v2_split"].eq(split)].copy().reset_index(drop=True)
    if result.empty:
        raise ValueError(f"Empty split: {split}")
    return result


def metrics_for(labels, predictions, probabilities) -> dict:
    labels = np.asarray(labels, dtype=int)
    predictions = np.asarray(predictions, dtype=int)
    probabilities = np.asarray(probabilities, dtype=float)
    result = {
        "accuracy": float(accuracy_score(labels, predictions)),
        "precision": float(precision_score(labels, predictions, zero_division=0)),
        "recall": float(recall_score(labels, predictions, zero_division=0)),
        "f1": float(f1_score(labels, predictions, zero_division=0)),
        "macro_f1": float(f1_score(labels, predictions, average="macro", zero_division=0)),
        "recall_class_0": float(recall_score(labels, predictions, labels=[0], average=None, zero_division=0)[0]),
        "recall_class_1": float(recall_score(labels, predictions, labels=[1], average=None, zero_division=0)[0]),
        "roc_auc": float(roc_auc_score(labels, probabilities)) if np.unique(labels).size == 2 else None,
        "pr_auc": float(average_precision_score(labels, probabilities)) if np.unique(labels).size == 2 else None,
        "confusion_matrix": confusion_matrix(labels, predictions, labels=[0, 1]).tolist(),
    }
    return result


class TextDataset(Dataset):
    def __init__(self, dataframe: pd.DataFrame, tokenizer):
        self.ids = dataframe["id"].astype(str).tolist()
        self.labels = torch.tensor(dataframe["label"].to_numpy(dtype=int), dtype=torch.long)
        self.encodings = tokenizer(
            dataframe["text"].fillna("").astype(str).tolist(),
            padding="max_length",
            truncation=True,
            max_length=MAX_LENGTH,
            return_tensors="pt",
        )

    def __len__(self):
        return len(self.labels)

    def __getitem__(self, index):
        item = {key: value[index] for key, value in self.encodings.items()}
        item["labels"] = self.labels[index]
        item["sample_index"] = torch.tensor(index, dtype=torch.long)
        return item


# END REGISTERED SOURCE BLOCK


In [99]:
%%project_source historical/v2/experiments/source_disjoint/run_source_disjoint.py 1
class ImageDataset(Dataset):
    def __init__(self, dataframe: pd.DataFrame, transform):
        self.df = dataframe.reset_index(drop=True)
        self.transform = transform

    def __len__(self):
        return len(self.df)

    def __getitem__(self, index):
        row = self.df.iloc[index]
        with Image.open(row["resolved_image_path"]) as image:
            tensor = self.transform(image.convert("RGB"))
        return {
            "image": tensor,
            "label": torch.tensor(int(row["label"]), dtype=torch.long),
            "sample_index": torch.tensor(index, dtype=torch.long),
        }


def image_transform():
    return transforms.Compose([
        transforms.Resize((224, 224)),
        transforms.ToTensor(),
        transforms.Normalize(mean=[0.485, 0.456, 0.406], std=[0.229, 0.224, 0.225]),
    ])


def worker_seed(worker_id: int) -> None:
    worker_seed_value = SEED + worker_id
    np.random.seed(worker_seed_value)
    random.seed(worker_seed_value)


def text_evaluate(model, loader, device):
    model.eval()
    labels, predictions, probabilities, indices = [], [], [], []
    total_loss = 0.0
    with torch.no_grad():
        for batch in loader:
            index = batch.pop("sample_index")
            cpu_labels = batch["labels"].numpy()
            batch = {key: value.to(device, non_blocking=True) for key, value in batch.items()}
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                output = model(**batch)
            probability = torch.softmax(output.logits, dim=1)[:, 1]
            prediction = (probability >= THRESHOLD).long()
            total_loss += float(output.loss.item())
            indices.extend(index.numpy().tolist())
            labels.extend(cpu_labels.tolist())
            predictions.extend(prediction.cpu().numpy().tolist())
            probabilities.extend(probability.cpu().float().numpy().tolist())
    result = metrics_for(labels, predictions, probabilities)
    result["loss"] = total_loss / len(loader)
    return result, np.asarray(indices), np.asarray(labels), np.asarray(predictions), np.asarray(probabilities)


def image_evaluate(model, loader, device):
    model.eval()
    labels, predictions, probabilities, indices = [], [], [], []
    total_loss = 0.0
    criterion = nn.CrossEntropyLoss()
    with torch.no_grad():
        for batch in loader:
            image = batch["image"].to(device, non_blocking=True)
            label = batch["label"].to(device, non_blocking=True)
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                logits = model(image)
                loss = criterion(logits, label)
            probability = torch.softmax(logits, dim=1)[:, 1]
            prediction = (probability >= THRESHOLD).long()
            total_loss += float(loss.item())
            indices.extend(batch["sample_index"].numpy().tolist())
            labels.extend(label.cpu().numpy().tolist())
            predictions.extend(prediction.cpu().numpy().tolist())
            probabilities.extend(probability.cpu().float().numpy().tolist())
    result = metrics_for(labels, predictions, probabilities)
    result["loss"] = total_loss / len(loader)
    return result, np.asarray(indices), np.asarray(labels), np.asarray(predictions), np.asarray(probabilities)


def prediction_frame(dataframe, indices, labels, predictions, probabilities, prefix: str) -> pd.DataFrame:
    indexed = dataframe.iloc[indices].reset_index(drop=True)
    if not np.array_equal(indexed["label"].to_numpy(dtype=int), labels):
        raise ValueError(f"Label alignment failed for {prefix}")
    return pd.DataFrame({
        "sample_id": indexed["id"].astype(str),
        "true_label": labels,
        f"{prefix}_probability_class1": probabilities,
        f"{prefix}_prediction": predictions,
    })


def stage_audit(root: Path) -> None:
    make_dirs(root)
    p = paths(root)
    if not SOURCE_MANIFEST.exists():
        raise FileNotFoundError(SOURCE_MANIFEST)
    if p["manifest"].exists():
        if hashlib.sha256(p["manifest"].read_bytes()).hexdigest() != hashlib.sha256(SOURCE_MANIFEST.read_bytes()).hexdigest():
            raise FileExistsError(f"An unrelated manifest already exists at {p['manifest']}")
    else:
        shutil.copy2(SOURCE_MANIFEST, p["manifest"])

    df = pd.read_parquet(p["manifest"])
    required = ["id", "label", "text", "image_path", "subreddit", "domain", "created_utc", "v2_split"]
    if list(df.columns) != required:
        raise ValueError(f"Unexpected schema: {df.columns.tolist()}")
    if df["id"].astype(str).duplicated().any():
        raise ValueError("Duplicate sample IDs")
    if set(df["v2_split"]) != {"train", "validation", "test"}:
        raise ValueError("Unexpected split labels")
    if set(df["label"].astype(int)) != {0, 1}:
        raise ValueError("Unexpected class labels")

    source_sets = {name: set(group["subreddit"].astype(str)) for name, group in df.groupby("v2_split")}
    overlap = {}
    names = sorted(source_sets)
    for i, left in enumerate(names):
        for right in names[i + 1:]:
            overlap[f"{left}__{right}"] = sorted(source_sets[left] & source_sets[right])
    if any(overlap.values()):
        raise ValueError(f"Source overlap found: {overlap}")

    records, unreadable, placeholders = [], [], []
    for row in df.itertuples(index=False):
        image_path = resolve_image_path(row.image_path)
        exists = image_path.is_file()
        readable = False
        digest = None
        error = None
        if exists:
            try:
                with Image.open(image_path) as image:
                    image.verify()
                readable = True
                digest = hashlib.sha256(image_path.read_bytes()).hexdigest()
            except Exception as exc:  # recorded in audit output
                error = repr(exc)
        if not readable:
            unreadable.append({"id": str(row.id), "path": str(image_path), "error": error or "missing"})
        if digest == PLACEHOLDER_SHA256:
            placeholders.append(str(row.id))
        records.append({"v2_split": row.v2_split, "label": int(row.label), "readable": readable})
    checks = pd.DataFrame(records)
    split_rows = []
    for split in ["train", "validation", "test"]:
        part = df[df["v2_split"].eq(split)]
        verified = checks[checks["v2_split"].eq(split)]
        split_rows.append({
            "split": split,
            "manifest_samples": int(len(part)),
            "retained_samples": int(verified["readable"].sum()),
            "removed_samples": int((~verified["readable"]).sum()),
            "removed_class_0": 0,
            "removed_class_1": 0,
            "class_0": int(part["label"].eq(0).sum()),
            "class_1": int(part["label"].eq(1).sum()),
            "class_1_rate": float(part["label"].mean()),
            "sources": int(part["subreddit"].nunique()),
        })
    if unreadable or placeholders:
        raise ValueError(f"Manifest contains {len(unreadable)} unreadable and {len(placeholders)} placeholder images")
    pd.DataFrame(split_rows).to_csv(p["manifests"] / "split_counts.csv", index=False)

    manifest_sha = hashlib.sha256(p["manifest"].read_bytes()).hexdigest()
    audit = {
        "source_manifest": str(SOURCE_MANIFEST),
        "isolated_manifest": str(p["manifest"]),
        "sha256": manifest_sha,
        "schema": {column: str(dtype) for column, dtype in df.dtypes.items()},
        "rows": int(len(df)),
        "duplicate_ids": 0,
        "blank_text": int(df["text"].fillna("").astype(str).str.strip().eq("").sum()),
        "source_overlap": overlap,
        "unreadable_images": unreadable,
        "known_placeholder_images": placeholders,
        "splits": split_rows,
        "positive_class": "1 (true)",
        "negative_class": "0 (fake or misleading)",
        "note": "The manifest was constructed from the existing cleaned multimodal pool, so its manifest and retained counts are equal.",
    }
    dump_json(p["audit"], audit)
    config = {
        "experiment": "source_disjoint",
        "created_utc": datetime.now(timezone.utc).isoformat(),
        "seed": SEED,
        "project_root": str(PROJECT_ROOT),
        "source_manifest": str(SOURCE_MANIFEST),
        "isolated_manifest": str(p["manifest"]),
        "manifest_sha256": manifest_sha,
        "split_counts": {row["split"]: row["retained_samples"] for row in split_rows},
        "positive_class": 1,
        "classification_threshold": THRESHOLD,
        "roberta": {"base_model": MODEL_NAME, "pretrained_base_weights": True, "max_length": MAX_LENGTH, "batch_size": 16, "optimizer": "AdamW", "learning_rate": 2e-5, "weight_decay": 0.01, "gradient_clipping": 1.0, "warmup_fraction": 0.10, "max_epochs": 3, "selection_metric": "validation_macro_f1", "checkpoint": str(p["roberta_checkpoint"])},
        "resnet50": {"base_model": "resnet50", "weights": "IMAGENET1K_V2", "fine_tune": "full network", "input_size": [224, 224], "batch_size": 32, "optimizer": "AdamW", "learning_rate": 1e-4, "weight_decay": 0.01, "max_epochs": 3, "selection_metric": "validation_macro_f1", "checkpoint": str(p["resnet_checkpoint"] / "best_model.pt")},
        "fusion": {"formula": "alpha * p_text + (1 - alpha) * p_image", "alpha_search": [round(x, 2) for x in np.arange(0, 1.0001, 0.05)], "selection_metric": "validation_macro_f1", "tie_break": "closest to 0.50, then lower alpha", "selected_alpha": None},
        "calibration": {"ece_bins": N_BINS, "convention": "confidence bins from 0.5 to 1.0"},
        "bootstrap": {"iterations": N_BOOTSTRAPS, "seed": SEED, "paired": True},
        "packages": {"python": platform.python_version(), "torch": torch.__version__, "torchvision": torchvision.__version__, "transformers": transformers.__version__, "pandas": pd.__version__, "numpy": np.__version__, "scikit_learn": sklearn.__version__, "scipy": scipy.__version__},
        "hardware": {"cuda_available": torch.cuda.is_available(), "cuda_version": torch.version.cuda, "gpu": torch.cuda.get_device_name(0) if torch.cuda.is_available() else None},
    }
    dump_json(p["config"], config)
    print(pd.DataFrame(split_rows).to_string(index=False))
    print(f"Audit saved: {p['audit']}")


# END REGISTERED SOURCE BLOCK


In [100]:
%%project_source historical/v2/experiments/source_disjoint/run_source_disjoint.py 2
def create_resnet() -> nn.Module:
    model = resnet50(weights=ResNet50_Weights.IMAGENET1K_V2)
    model.fc = nn.Linear(model.fc.in_features, 2)
    return model


def stage_smoke(root: Path) -> None:
    set_seed()
    df = load_manifest(root)
    train = split_df(df, "train").sample(n=32, random_state=SEED).reset_index(drop=True)
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    tokenizer = AutoTokenizer.from_pretrained(MODEL_NAME)
    text_loader = DataLoader(TextDataset(train, tokenizer), batch_size=8, shuffle=False)
    text_model = AutoModelForSequenceClassification.from_pretrained(MODEL_NAME, num_labels=2).to(device)
    text_batch = next(iter(text_loader))
    text_indices = text_batch.pop("sample_index")
    with torch.no_grad(), torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
        text_out = text_model(**{key: value.to(device) for key, value in text_batch.items()})
    image_loader = DataLoader(ImageDataset(train, image_transform()), batch_size=4, shuffle=False, num_workers=0)
    image_model = create_resnet().to(device)
    image_batch = next(iter(image_loader))
    with torch.no_grad(), torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
        image_logits = image_model(image_batch["image"].to(device))
    if text_out.logits.shape != (8, 2) or image_logits.shape != (4, 2):
        raise ValueError("Unexpected smoke-test output shape")
    if not np.array_equal(text_batch["labels"].numpy(), train.iloc[text_indices.numpy()]["label"].to_numpy()):
        raise ValueError("Text labels are not aligned")
    if not np.array_equal(image_batch["label"].numpy(), train.iloc[image_batch["sample_index"].numpy()]["label"].to_numpy()):
        raise ValueError("Image labels are not aligned")
    result = {"passed": True, "device": str(device), "gpu": torch.cuda.get_device_name(0) if device.type == "cuda" else None, "text_batch_shape": list(text_out.logits.shape), "image_batch_shape": list(image_logits.shape), "labels_aligned": True, "output_root": str(root)}
    dump_json(paths(root)["logs"] / "smoke_test.json", result)
    print(json.dumps(result, indent=2))


def train_roberta(root: Path, epochs: int, batch_size: int) -> None:
    p = paths(root)
    if (p["roberta_checkpoint"] / "model.safetensors").exists() or (p["roberta_checkpoint"] / "pytorch_model.bin").exists():
        raise FileExistsError("RoBERTa checkpoint already exists; refusing to overwrite it")
    set_seed()
    df = load_manifest(root)
    train, validation = split_df(df, "train"), split_df(df, "validation")
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    tokenizer = AutoTokenizer.from_pretrained(MODEL_NAME)
    train_loader = DataLoader(TextDataset(train, tokenizer), batch_size=batch_size, shuffle=True, num_workers=0, pin_memory=device.type == "cuda", generator=torch.Generator().manual_seed(SEED))
    validation_loader = DataLoader(TextDataset(validation, tokenizer), batch_size=batch_size, shuffle=False, num_workers=0, pin_memory=device.type == "cuda")
    model = AutoModelForSequenceClassification.from_pretrained(MODEL_NAME, num_labels=2).to(device)
    optimizer = AdamW(model.parameters(), lr=2e-5, weight_decay=0.01)
    total_steps = len(train_loader) * epochs
    scheduler = get_linear_schedule_with_warmup(optimizer, num_warmup_steps=int(total_steps * 0.10), num_training_steps=total_steps)
    scaler = torch.amp.GradScaler("cuda", enabled=device.type == "cuda")
    history, best = [], -1.0
    for epoch in range(1, epochs + 1):
        model.train()
        total_loss = 0.0
        for step, batch in enumerate(train_loader, 1):
            batch.pop("sample_index")
            batch = {key: value.to(device, non_blocking=True) for key, value in batch.items()}
            optimizer.zero_grad(set_to_none=True)
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                output = model(**batch)
                loss = output.loss
            scaler.scale(loss).backward()
            scaler.unscale_(optimizer)
            torch.nn.utils.clip_grad_norm_(model.parameters(), 1.0)
            scaler.step(optimizer)
            scaler.update()
            scheduler.step()
            total_loss += float(loss.item())
            if step % 100 == 0:
                print(f"RoBERTa epoch {epoch} step {step}/{len(train_loader)} loss={total_loss/step:.4f}", flush=True)
        val_metrics, indices, labels, preds, probs = text_evaluate(model, validation_loader, device)
        record = {"epoch": epoch, "train_loss": total_loss / len(train_loader), **{f"validation_{k}": v for k, v in val_metrics.items() if k != "confusion_matrix"}}
        history.append(record)
        print(json.dumps(record, allow_nan=False), flush=True)
        if val_metrics["macro_f1"] > best:
            best = val_metrics["macro_f1"]
            model.save_pretrained(p["roberta_checkpoint"])
            tokenizer.save_pretrained(p["roberta_checkpoint"])
            prediction_frame(validation, indices, labels, preds, probs, "roberta").to_csv(p["predictions"] / "roberta_validation.csv", index=False)
            dump_json(p["metrics"] / "roberta_best_validation.json", {"best_epoch": epoch, "metrics": val_metrics, "checkpoint": str(p["roberta_checkpoint"])})
    pd.DataFrame(history).to_csv(p["metrics"] / "roberta_training_history.csv", index=False)
    print(f"Best validation macro F1: {best:.6f}")


def train_resnet(root: Path, epochs: int, batch_size: int, num_workers: int) -> None:
    p = paths(root)
    checkpoint_path = p["resnet_checkpoint"] / "best_model.pt"
    if checkpoint_path.exists():
        raise FileExistsError("ResNet checkpoint already exists; refusing to overwrite it")
    set_seed()
    df = load_manifest(root)
    train, validation = split_df(df, "train"), split_df(df, "validation")
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")
    loader_args = {"num_workers": num_workers, "pin_memory": device.type == "cuda", "worker_init_fn": worker_seed}
    if num_workers > 0:
        loader_args["persistent_workers"] = True
    train_loader = DataLoader(ImageDataset(train, image_transform()), batch_size=batch_size, shuffle=True, generator=torch.Generator().manual_seed(SEED), **loader_args)
    validation_loader = DataLoader(ImageDataset(validation, image_transform()), batch_size=batch_size, shuffle=False, **loader_args)
    model = create_resnet().to(device)
    criterion = nn.CrossEntropyLoss()
    optimizer = AdamW(model.parameters(), lr=1e-4, weight_decay=0.01)
    scaler = torch.amp.GradScaler("cuda", enabled=device.type == "cuda")
    history, best = [], -1.0
    for epoch in range(1, epochs + 1):
        model.train()
        total_loss = 0.0
        for step, batch in enumerate(train_loader, 1):
            images = batch["image"].to(device, non_blocking=True)
            labels = batch["label"].to(device, non_blocking=True)
            optimizer.zero_grad(set_to_none=True)
            with torch.autocast(device_type="cuda", dtype=torch.float16, enabled=device.type == "cuda"):
                logits = model(images)
                loss = criterion(logits, labels)
            scaler.scale(loss).backward()
            scaler.unscale_(optimizer)
            torch.nn.utils.clip_grad_norm_(model.parameters(), 1.0)
            scaler.step(optimizer)
            scaler.update()
            total_loss += float(loss.item())
            if step % 50 == 0:
                print(f"ResNet epoch {epoch} step {step}/{len(train_loader)} loss={total_loss/step:.4f}", flush=True)
        val_metrics, indices, labels, preds, probs = image_evaluate(model, validation_loader, device)
        record = {"epoch": epoch, "train_loss": total_loss / len(train_loader), **{f"validation_{k}": v for k, v in val_metrics.items() if k != "confusion_matrix"}}
        history.append(record)
        print(json.dumps(record, allow_nan=False), flush=True)
        if val_metrics["macro_f1"] > best:
            best = val_metrics["macro_f1"]
            torch.save({"model_state_dict": model.state_dict(), "model": "resnet50", "weights": "IMAGENET1K_V2", "num_classes": 2, "best_epoch": epoch, "validation_macro_f1": best}, checkpoint_path)
            prediction_frame(validation, indices, labels, preds, probs, "resnet").to_csv(p["predictions"] / "resnet_validation.csv", index=False)
            dump_json(p["metrics"] / "resnet_best_validation.json", {"best_epoch": epoch, "metrics": val_metrics, "checkpoint": str(checkpoint_path)})
    pd.DataFrame(history).to_csv(p["metrics"] / "resnet_training_history.csv", index=False)
    print(f"Best validation macro F1: {best:.6f}")


def stage_lock(root: Path) -> None:
    p = paths(root)
    if p["lock"].exists():
        raise FileExistsError("Validation lock already exists; refusing to replace it")
    text = pd.read_csv(p["predictions"] / "roberta_validation.csv")
    image = pd.read_csv(p["predictions"] / "resnet_validation.csv")
    merged = text.merge(image, on=["sample_id", "true_label"], validate="one_to_one")
    expected = len(split_df(load_manifest(root), "validation"))
    if len(merged) != expected:
        raise ValueError(f"Paired validation count {len(merged)} does not equal {expected}")
    merged.to_csv(p["predictions"] / "validation_predictions.csv", index=False)
    rows = []
    y = merged["true_label"].to_numpy(dtype=int)
    for alpha in np.arange(0, 1.0001, 0.05):
        probability = alpha * merged["roberta_probability_class1"].to_numpy() + (1 - alpha) * merged["resnet_probability_class1"].to_numpy()
        pred = (probability >= THRESHOLD).astype(int)
        score = metrics_for(y, pred, probability)
        rows.append({"alpha_text": round(float(alpha), 2), "alpha_image": round(float(1-alpha), 2), **{k: v for k, v in score.items() if k not in {"confusion_matrix", "recall_class_0", "recall_class_1"}}})
    search = pd.DataFrame(rows)
    search.to_csv(p["metrics"] / "validation_alpha_search.csv", index=False)
    maximum = search["macro_f1"].max()
    tied = search[np.isclose(search["macro_f1"], maximum)].copy()
    tied["distance_from_half"] = (tied["alpha_text"] - 0.5).abs()
    selected = tied.sort_values(["distance_from_half", "alpha_text"], ascending=[True, True]).iloc[0]

    # Optional fair text control: tune threshold and Platt calibration on validation only.
    threshold_rows = []
    for threshold in np.arange(0.05, 0.951, 0.01):
        pred = (merged["roberta_probability_class1"].to_numpy() >= threshold).astype(int)
        threshold_rows.append({"threshold": round(float(threshold), 2), "macro_f1": f1_score(y, pred, average="macro", zero_division=0)})
    threshold_search = pd.DataFrame(threshold_rows)
    threshold_search.to_csv(p["metrics"] / "roberta_validation_threshold_search.csv", index=False)
    threshold_best = threshold_search.sort_values(["macro_f1", "threshold"], ascending=[False, True]).iloc[0]
    calibrator = LogisticRegression(random_state=SEED).fit(merged[["roberta_probability_class1"]], y)
    dump_json(p["metrics"] / "fair_text_validation_control.json", {"selected_threshold": float(threshold_best["threshold"]), "validation_macro_f1": float(threshold_best["macro_f1"]), "platt_coefficient": float(calibrator.coef_[0, 0]), "platt_intercept": float(calibrator.intercept_[0])})

    lock = {"locked_utc": datetime.now(timezone.utc).isoformat(), "selection_partition": "validation", "paired_validation_samples": int(len(merged)), "selection_metric": "macro_f1", "selected_alpha_text": float(selected["alpha_text"]), "selected_alpha_image": float(selected["alpha_image"]), "validation_macro_f1": float(selected["macro_f1"]), "classification_threshold": THRESHOLD, "tied_alpha_values": tied["alpha_text"].astype(float).tolist(), "tie_break": "closest to 0.50, then lower alpha", "roberta_checkpoint": str(p["roberta_checkpoint"]), "resnet_checkpoint": str(p["resnet_checkpoint"] / "best_model.pt")}
    dump_json(p["lock"], lock)
    config = json.loads(p["config"].read_text(encoding="utf-8"))
    config["fusion"]["selected_alpha"] = lock["selected_alpha_text"]
    config["fusion"]["locked_utc"] = lock["locked_utc"]
    dump_json(p["config"], config)
    print(json.dumps(lock, indent=2))


# END REGISTERED SOURCE BLOCK


In [101]:
%%project_source historical/v2/experiments/source_disjoint/run_source_disjoint.py 3
def ece(labels, probabilities, n_bins=N_BINS):
    labels = np.asarray(labels, dtype=int)
    probabilities = np.asarray(probabilities, dtype=float)
    predictions = (probabilities >= 0.5).astype(int)
    confidence = np.maximum(probabilities, 1 - probabilities)
    correctness = (predictions == labels).astype(float)
    edges = np.linspace(0.5, 1.0, n_bins + 1)
    value, rows = 0.0, []
    for index, (lower, upper) in enumerate(zip(edges[:-1], edges[1:])):
        mask = (confidence >= lower) & (confidence <= upper if index == n_bins - 1 else confidence < upper)
        count = int(mask.sum())
        mean_confidence = float(confidence[mask].mean()) if count else None
        accuracy = float(correctness[mask].mean()) if count else None
        gap = abs(accuracy - mean_confidence) if count else None
        if count:
            value += count / len(labels) * gap
        rows.append({"bin_lower": float(lower), "bin_upper": float(upper), "count": count, "mean_confidence": mean_confidence, "accuracy": accuracy, "gap": gap})
    return float(value), rows


def calibration_for(name, labels, probabilities):
    clipped = np.clip(np.asarray(probabilities, dtype=float), 1e-7, 1 - 1e-7)
    ece_value, bins = ece(labels, clipped)
    return {"model": name, "brier": float(brier_score_loss(labels, clipped)), "log_loss": float(log_loss(labels, clipped)), "ece": ece_value}, bins


def bootstrap(root: Path, y, models: dict[str, tuple[np.ndarray, np.ndarray]]) -> pd.DataFrame:
    rng = np.random.default_rng(SEED)
    text_pred, text_prob = models["roberta"]
    fusion_pred, fusion_prob = models["late_fusion"]
    observed_text = metrics_for(y, text_pred, text_prob)
    observed_fusion = metrics_for(y, fusion_pred, fusion_prob)
    names = ["accuracy", "f1", "macro_f1", "roc_auc", "pr_auc"]
    values = {name: [] for name in names}
    for _ in range(N_BOOTSTRAPS):
        idx = rng.integers(0, len(y), size=len(y))
        ys = y[idx]
        basic_text = metrics_for(ys, text_pred[idx], text_prob[idx])
        basic_fusion = metrics_for(ys, fusion_pred[idx], fusion_prob[idx])
        for name in names:
            if basic_text[name] is not None and basic_fusion[name] is not None:
                values[name].append(basic_fusion[name] - basic_text[name])
    pd.DataFrame({name: pd.Series(series) for name, series in values.items()}).to_csv(paths(root)["bootstrap"] / "paired_differences.csv", index=False)
    rows = []
    for name in names:
        series = np.asarray(values[name])
        rows.append({"metric": name, "difference": observed_fusion[name] - observed_text[name], "ci_lower": float(np.percentile(series, 2.5)), "ci_upper": float(np.percentile(series, 97.5)), "valid_iterations": int(len(series)), "requested_iterations": N_BOOTSTRAPS})
    result = pd.DataFrame(rows)
    result.to_csv(paths(root)["metrics"] / "statistical_comparison.csv", index=False)
    return result


def reliability_plot(root: Path, bins_by_model: dict[str, list[dict]]) -> None:
    fig, ax = plt.subplots(figsize=(7, 6))
    ax.plot([0.5, 1.0], [0.5, 1.0], color="black", linestyle=":", label="Perfect calibration")
    for name, rows in bins_by_model.items():
        frame = pd.DataFrame(rows).dropna(subset=["mean_confidence", "accuracy"])
        ax.plot(frame["mean_confidence"], frame["accuracy"], marker="o", label=name)
    ax.set(xlabel="Mean confidence", ylabel="Observed accuracy", xlim=(0.5, 1.0), ylim=(0.5, 1.0), title="Source-disjoint test reliability")
    ax.legend()
    fig.tight_layout()
    fig.savefig(paths(root)["figures"] / "reliability_diagram.png", dpi=180)
    plt.close(fig)


def markdown_table(frame: pd.DataFrame, decimals: int = 4) -> str:
    """Render a small DataFrame without the optional tabulate dependency."""
    display = frame.copy()
    for column in display.select_dtypes(include=["float", "floating"]).columns:
        display[column] = display[column].map(lambda value: "" if pd.isna(value) else f"{value:.{decimals}f}")
    headers = [str(column) for column in display.columns]
    lines = ["| " + " | ".join(headers) + " |", "| " + " | ".join(["---"] * len(headers)) + " |"]
    for row in display.itertuples(index=False, name=None):
        lines.append("| " + " | ".join(str(value).replace("|", "\\|") for value in row) + " |")
    return "\n".join(lines)


def stage_test(root: Path, text_batch: int, image_batch: int, num_workers: int) -> None:
    p = paths(root)
    final_predictions_path = p["predictions"] / "test_predictions.csv"
    if final_predictions_path.exists():
        raise FileExistsError("Test predictions already exist; refusing to evaluate the locked test twice")
    lock = json.loads(p["lock"].read_text(encoding="utf-8"))
    alpha = float(lock["selected_alpha_text"])
    set_seed()
    test = split_df(load_manifest(root), "test")
    device = torch.device("cuda" if torch.cuda.is_available() else "cpu")

    tokenizer = AutoTokenizer.from_pretrained(p["roberta_checkpoint"])
    text_loader = DataLoader(TextDataset(test, tokenizer), batch_size=text_batch, shuffle=False, num_workers=0, pin_memory=device.type == "cuda")
    text_model = AutoModelForSequenceClassification.from_pretrained(p["roberta_checkpoint"]).to(device)
    _, ti, ty, tp, tprob = text_evaluate(text_model, text_loader, device)
    text_frame = prediction_frame(test, ti, ty, tp, tprob, "roberta")
    del text_model
    if device.type == "cuda":
        torch.cuda.empty_cache()

    loader_args = {"num_workers": num_workers, "pin_memory": device.type == "cuda", "worker_init_fn": worker_seed}
    if num_workers > 0:
        loader_args["persistent_workers"] = True
    image_loader = DataLoader(ImageDataset(test, image_transform()), batch_size=image_batch, shuffle=False, **loader_args)
    image_model = create_resnet().to(device)
    checkpoint = torch.load(p["resnet_checkpoint"] / "best_model.pt", map_location=device, weights_only=True)
    image_model.load_state_dict(checkpoint["model_state_dict"])
    _, ii, iy, ip, iprob = image_evaluate(image_model, image_loader, device)
    image_frame = prediction_frame(test, ii, iy, ip, iprob, "resnet")

    predictions = text_frame.merge(image_frame, on=["sample_id", "true_label"], validate="one_to_one")
    diagnostics = test[["id", "subreddit"]].rename(columns={"id": "sample_id"})
    predictions = predictions.merge(diagnostics, on="sample_id", validate="one_to_one")
    predictions["fusion_probability_class1"] = alpha * predictions["roberta_probability_class1"] + (1 - alpha) * predictions["resnet_probability_class1"]
    predictions["fusion_prediction"] = (predictions["fusion_probability_class1"] >= THRESHOLD).astype(int)
    predictions.to_csv(final_predictions_path, index=False)

    y = predictions["true_label"].to_numpy(dtype=int)
    model_arrays = {
        "roberta": (predictions["roberta_prediction"].to_numpy(dtype=int), predictions["roberta_probability_class1"].to_numpy()),
        "resnet50": (predictions["resnet_prediction"].to_numpy(dtype=int), predictions["resnet_probability_class1"].to_numpy()),
        "late_fusion": (predictions["fusion_prediction"].to_numpy(dtype=int), predictions["fusion_probability_class1"].to_numpy()),
    }
    metric_rows, full_metrics = [], {}
    calibration_rows, bins_by_model = [], {}
    for name, (pred, prob) in model_arrays.items():
        values = metrics_for(y, pred, prob)
        full_metrics[name] = values
        cal, bins = calibration_for(name, y, prob)
        calibration_rows.append(cal)
        bins_by_model[name] = bins
        pd.DataFrame(bins).to_csv(p["calibration"] / f"{name}_bins.csv", index=False)
        metric_rows.append({"model": name, **{key: value for key, value in values.items() if key != "confusion_matrix"}, **{key: value for key, value in cal.items() if key != "model"}})
    metric_summary = pd.DataFrame(metric_rows)
    metric_summary.to_csv(p["metrics"] / "summary.csv", index=False)
    dump_json(p["metrics"] / "summary.json", {"test_samples": len(predictions), "selected_alpha_text": alpha, "models": full_metrics})
    calibration_frame = pd.DataFrame(calibration_rows)
    calibration_frame.to_csv(p["calibration"] / "calibration_metrics.csv", index=False)
    dump_json(p["calibration"] / "calibration_metrics.json", {"n_bins": N_BINS, "convention": "confidence bins from 0.5 to 1.0", "models": calibration_rows})
    reliability_plot(root, bins_by_model)

    cr = model_arrays["roberta"][0] == y
    ci = model_arrays["resnet50"][0] == y
    cf = model_arrays["late_fusion"][0] == y
    b = int(np.sum(cr & ~cf))
    c = int(np.sum(~cr & cf))
    mcnemar_p = float(binomtest(min(b, c), n=b + c, p=0.5, alternative="two-sided").pvalue) if b + c else 1.0
    mcnemar = {"both_correct": int(np.sum(cr & cf)), "both_wrong": int(np.sum(~cr & ~cf)), "roberta_correct_fusion_wrong": b, "fusion_correct_roberta_wrong": c, "discordant": b + c, "exact_p_value": mcnemar_p}
    dump_json(p["metrics"] / "mcnemar.json", mcnemar)
    stats = bootstrap(root, y, model_arrays)
    complementarity = {
        "roberta_vs_fusion": mcnemar,
        "roberta_vs_resnet_disagreements": int(np.sum(model_arrays["roberta"][0] != model_arrays["resnet50"][0])),
        "roberta_only_correct": int(np.sum(cr & ~ci)),
        "resnet_only_correct": int(np.sum(~cr & ci)),
        "image_correct_text_wrong_recovered_by_fusion": int(np.sum(~cr & ci & cf)),
        "text_correct_image_wrong_preserved_by_fusion": int(np.sum(cr & ~ci & cf)),
    }
    dump_json(p["metrics"] / "error_complementarity.json", complementarity)

    # Apply the validation-selected fair text threshold and Platt model once to test.
    fair = json.loads((p["metrics"] / "fair_text_validation_control.json").read_text(encoding="utf-8"))
    tuned_pred = (model_arrays["roberta"][1] >= fair["selected_threshold"]).astype(int)
    z = fair["platt_intercept"] + fair["platt_coefficient"] * model_arrays["roberta"][1]
    platt_prob = 1 / (1 + np.exp(-z))
    pd.DataFrame([
        {"control": "validation_tuned_threshold", "threshold": fair["selected_threshold"], **{k: v for k, v in metrics_for(y, tuned_pred, model_arrays["roberta"][1]).items() if k != "confusion_matrix"}},
        {"control": "validation_platt_calibration", "threshold": 0.5, **{k: v for k, v in metrics_for(y, (platt_prob >= 0.5).astype(int), platt_prob).items() if k != "confusion_matrix"}},
    ]).to_csv(p["metrics"] / "fair_text_test_control.csv", index=False)

    original = {"roberta": {"accuracy": 0.8046, "macro_f1": 0.8000, "roc_auc": 0.8846, "pr_auc": 0.9027}, "resnet50": {"accuracy": 0.7382, "macro_f1": 0.7275, "roc_auc": 0.7976, "pr_auc": 0.8053}, "late_fusion": {"accuracy": 0.8242, "macro_f1": 0.8188, "roc_auc": 0.8993, "pr_auc": 0.9097}}
    penalty_rows = []
    for name in original:
        for metric, old in original[name].items():
            penalty_rows.append({"model": name, "metric": metric, "ordinary_locked_holdout": old, "source_disjoint": full_metrics[name][metric], "change_source_disjoint_minus_ordinary": full_metrics[name][metric] - old})
    pd.DataFrame(penalty_rows).to_csv(p["metrics"] / "generalisation_penalty.csv", index=False)

    counts = pd.read_csv(p["manifests"] / "split_counts.csv")
    macro_row = stats[stats["metric"].eq("macro_f1")].iloc[0]
    best_text = json.loads((p["metrics"] / "roberta_best_validation.json").read_text(encoding="utf-8"))
    best_image = json.loads((p["metrics"] / "resnet_best_validation.json").read_text(encoding="utf-8"))
    lines = [
        "# Source-disjoint evaluation results", "",
        "## Dataset and split verification", "",
        "The manifest assigns every subreddit to one partition. No subreddit appears in more than one split. Both labels occur in every split. All image files opened correctly and the known regional-unavailable placeholder was absent.", "",
        markdown_table(counts), "",
        "The source-disjoint manifest was created from the existing cleaned multimodal pool. The manifest count is therefore also the final usable count, with no further removals in this run.", "",
        "## Locked validation choices", "",
        f"RoBERTa checkpoint: `{best_text['checkpoint']}` (epoch {best_text['best_epoch']}).", "",
        f"ResNet-50 checkpoint: `{best_image['checkpoint']}` (epoch {best_image['best_epoch']}).", "",
        f"Validation selected alpha = {alpha:.2f} for RoBERTa and {1-alpha:.2f} for ResNet-50. The classification threshold remained 0.50.", "",
        "The complete search is in `metrics/validation_alpha_search.csv`.", "",
        "## Source-disjoint test performance", "", markdown_table(metric_summary), "",
        "## Calibration", "", markdown_table(calibration_frame), "",
        "Lower Brier score, log loss and ECE indicate better calibration.", "",
        "## Paired statistical comparison", "",
        f"Late fusion and RoBERTa were compared on {len(y):,} paired test cases. Both were correct on {mcnemar['both_correct']:,}; both were wrong on {mcnemar['both_wrong']:,}. RoBERTa alone was correct on {b:,} and fusion alone on {c:,}. The exact McNemar p-value was {mcnemar_p:.6g}.", "",
        markdown_table(stats), "",
        "## Error complementarity", "",
        f"RoBERTa and ResNet-50 disagreed on {complementarity['roberta_vs_resnet_disagreements']:,} cases. RoBERTa alone was correct on {complementarity['roberta_only_correct']:,}; ResNet-50 alone was correct on {complementarity['resnet_only_correct']:,}. Late fusion recovered {complementarity['image_correct_text_wrong_recovered_by_fusion']:,} image-correct/text-wrong cases and preserved {complementarity['text_correct_image_wrong_preserved_by_fusion']:,} text-correct/image-wrong cases.", "",
        "## Interpretation", "",
        f"Removing subreddit overlap changed RoBERTa macro F1 by {full_metrics['roberta']['macro_f1']-0.8000:+.4f}, ResNet-50 by {full_metrics['resnet50']['macro_f1']-0.7275:+.4f}, and late fusion by {full_metrics['late_fusion']['macro_f1']-0.8188:+.4f} compared with the ordinary locked holdout. Late fusion changed macro F1 over RoBERTa by {full_metrics['late_fusion']['macro_f1']-full_metrics['roberta']['macro_f1']:+.4f}. Its paired 95% bootstrap interval was [{macro_row['ci_lower']:+.4f}, {macro_row['ci_upper']:+.4f}]. Validation selected zero text weight, so the locked late-fusion result is identical to ResNet-50 and does not show a benefit from combining modalities. These figures measure transfer to unseen subreddit groups rather than performance on the earlier mixed-source holdout.", "",
    ]
    (p["reports"] / "source_disjoint_results.md").write_text("\n".join(lines), encoding="utf-8")
    config = json.loads(p["config"].read_text(encoding="utf-8"))
    config["test_evaluated_utc"] = datetime.now(timezone.utc).isoformat()
    config["test_predictions"] = str(final_predictions_path)
    dump_json(p["config"], config)
    print(metric_summary.to_string(index=False))
    print(json.dumps(mcnemar, indent=2))


# END REGISTERED SOURCE BLOCK


In [102]:
%%project_source historical/v2/experiments/source_disjoint/run_source_disjoint.py 4
def main() -> None:
    parser = argparse.ArgumentParser()
    parser.add_argument("stage", choices=["audit", "smoke", "train-roberta", "train-resnet", "lock", "test"])
    parser.add_argument("--experiment-root", type=Path, default=DEFAULT_EXPERIMENT_ROOT)
    parser.add_argument("--epochs", type=int, default=3)
    parser.add_argument("--batch-size", type=int)
    parser.add_argument("--num-workers", type=int, default=2)
    args = parser.parse_args()
    root = args.experiment_root.resolve()
    if args.stage == "audit": stage_audit(root)
    elif args.stage == "smoke": stage_smoke(root)
    elif args.stage == "train-roberta": train_roberta(root, args.epochs, args.batch_size or 16)
    elif args.stage == "train-resnet": train_resnet(root, args.epochs, args.batch_size or 32, args.num_workers)
    elif args.stage == "lock": stage_lock(root)
    elif args.stage == "test": stage_test(root, args.batch_size or 16, 32, args.num_workers)


if __name__ == "__main__":
    main()
# END REGISTERED SOURCE BLOCK


#### Earlier local file: `v2/experiments/source_disjoint/build_report.py`

In [103]:
%%project_source historical/v2/experiments/source_disjoint/build_report.py 0
"""Build the source-disjoint Markdown report from already saved outputs."""
from __future__ import annotations

import json
from datetime import datetime, timezone
from pathlib import Path

import pandas as pd


ROOT = Path(r"F:\data sci\project\v2\experiments\source_disjoint")


def table(frame: pd.DataFrame, decimals: int = 4) -> str:
    data = frame.copy()
    for column in data.select_dtypes(include=["float", "floating"]).columns:
        data[column] = data[column].map(lambda value: "" if pd.isna(value) else f"{value:.{decimals}f}")
    lines = [
        "| " + " | ".join(map(str, data.columns)) + " |",
        "| " + " | ".join(["---"] * len(data.columns)) + " |",
    ]
    for row in data.itertuples(index=False, name=None):
        lines.append("| " + " | ".join(str(value).replace("|", "\\|") for value in row) + " |")
    return "\n".join(lines)


def load_json(relative: str):
    return json.loads((ROOT / relative).read_text(encoding="utf-8"))


counts = pd.read_csv(ROOT / "manifests/split_counts.csv")
summary = pd.read_csv(ROOT / "metrics/summary.csv")
calibration = pd.read_csv(ROOT / "calibration/calibration_metrics.csv")
stats = pd.read_csv(ROOT / "metrics/statistical_comparison.csv")
alpha_search = pd.read_csv(ROOT / "metrics/validation_alpha_search.csv")
penalty = pd.read_csv(ROOT / "metrics/generalisation_penalty.csv")
lock = load_json("metrics/validation_lock.json")
mcnemar = load_json("metrics/mcnemar.json")
errors = load_json("metrics/error_complementarity.json")
text_best = load_json("metrics/roberta_best_validation.json")
image_best = load_json("metrics/resnet_best_validation.json")

metrics = summary.set_index("model")
macro = stats.set_index("metric").loc["macro_f1"]
alpha = lock["selected_alpha_text"]

lines = [
    "# Source-disjoint evaluation results",
    "",
    "## Dataset and split verification",
    "",
    "The copied manifest contains 17,056 cleaned multimodal samples. Each subreddit belongs to one partition only and both labels appear in each split. All image paths resolve, every image opens correctly and the regional-unavailable placeholder is absent. Sample IDs are unique and all text fields are non-empty.",
    "",
    table(counts),
    "",
    "The source-disjoint manifest was built from the existing cleaned multimodal pool. Its manifest count is also its final usable count, so this run removed no further samples from either class.",
    "",
    "## Training and locked validation choices",
    "",
    "RoBERTa-base and ResNet-50 were trained from their pretrained base weights using only the source-disjoint training split. Subreddit, domain, timestamp and engagement fields were not model inputs. Both models used a maximum of three epochs and the best checkpoint was chosen by validation macro F1.",
    "",
    f"RoBERTa checkpoint: `{text_best['checkpoint']}`. Epoch {text_best['best_epoch']} was selected with validation macro F1 {text_best['metrics']['macro_f1']:.4f}.",
    "",
    f"ResNet-50 checkpoint: `{image_best['checkpoint']}`. Epoch {image_best['best_epoch']} was selected with validation macro F1 {image_best['metrics']['macro_f1']:.4f}.",
    "",
    f"The validation search selected α = {alpha:.2f} for RoBERTa and {1-alpha:.2f} for ResNet-50 at threshold 0.50. There was no tie. Since α is zero, the locked late-fusion model is numerically identical to ResNet-50. It should not be described as a benefit from combining modalities.",
    "",
    "The full 21-point search is saved in `metrics/validation_alpha_search.csv`.",
    "",
    "## Source-disjoint test performance",
    "",
    table(summary),
    "",
    "RoBERTa remained the stronger unimodal model on the three unseen test subreddits. ResNet-50 retained predictive information but scored below RoBERTa. The validation-selected late fusion also scored below RoBERTa because validation assigned zero weight to text.",
    "",
    "## Calibration",
    "",
    table(calibration),
    "",
    "ResNet-50 and the locked fusion had lower ECE, while RoBERTa had lower Brier score and log loss. ECE uses the project convention of ten confidence bins from 0.5 to 1.0.",
    "",
    "## McNemar test",
    "",
    f"Both RoBERTa and fusion were correct on {mcnemar['both_correct']:,} cases and both were wrong on {mcnemar['both_wrong']:,}. RoBERTa alone was correct on {mcnemar['roberta_correct_fusion_wrong']:,}; fusion alone was correct on {mcnemar['fusion_correct_roberta_wrong']:,}. The exact two-sided McNemar p-value was {mcnemar['exact_p_value']:.6g}.",
    "",
    "The direction favours RoBERTa because it won more discordant cases.",
    "",
    "## Paired bootstrap confidence intervals",
    "",
    table(stats),
    "",
    f"The fusion-minus-RoBERTa macro F1 difference was {macro['difference']:+.4f}, with a 95% paired bootstrap interval of [{macro['ci_lower']:+.4f}, {macro['ci_upper']:+.4f}]. The interval does not cross zero and favours RoBERTa.",
    "",
    "## Error complementarity",
    "",
    f"RoBERTa and ResNet-50 disagreed on {errors['roberta_vs_resnet_disagreements']:,} test cases. RoBERTa alone was correct on {errors['roberta_only_correct']:,}; ResNet-50 alone was correct on {errors['resnet_only_correct']:,}. The locked fusion recovered all {errors['image_correct_text_wrong_recovered_by_fusion']:,} image-correct/text-wrong cases because it equals the image model, but it preserved none of the {errors['roberta_only_correct']:,} text-correct/image-wrong cases.",
    "",
    "The disagreement count shows that the modalities make different errors. The selected coefficient did not use that complementarity on test because the two validation subreddits favoured an image-only decision.",
    "",
    "## Change from the ordinary locked holdout",
    "",
    table(penalty),
    "",
    f"RoBERTa macro F1 fell from 0.8000 to {metrics.loc['roberta', 'macro_f1']:.4f}, a change of {metrics.loc['roberta', 'macro_f1']-0.8000:+.4f}. ResNet-50 fell from 0.7275 to {metrics.loc['resnet50', 'macro_f1']:.4f}, a change of {metrics.loc['resnet50', 'macro_f1']-0.7275:+.4f}. Locked late fusion fell from 0.8188 to {metrics.loc['late_fusion', 'macro_f1']:.4f}, a change of {metrics.loc['late_fusion', 'macro_f1']-0.8188:+.4f}.",
    "",
    "## Interpretation",
    "",
    "Removing source overlap produced a clear generalisation penalty for all three reported systems. RoBERTa still transferred better than ResNet-50 on the test sources. The image model retained useful signal, shown by its ROC AUC and the cases it alone classified correctly.",
    "",
    "Late fusion did not outperform RoBERTa in this experiment. Its validation-selected coefficient removed the text contribution, then underperformed RoBERTa on test by 0.0825 macro F1. The confidence interval and McNemar result support that direction. This also exposes a limit in the split: validation contains only two subreddits and test contains three. Model and fusion selection can depend heavily on which whole sources enter each partition. The result is still useful because it shows how performance and modality weighting change when source overlap is removed.",
    "",
]

report_path = ROOT / "reports/source_disjoint_results.md"
report_path.parent.mkdir(parents=True, exist_ok=True)
report_path.write_text("\n".join(lines), encoding="utf-8")

config_path = ROOT / "experiment_config.json"
config = json.loads(config_path.read_text(encoding="utf-8"))
config["test_evaluated_utc"] = datetime.now(timezone.utc).isoformat()
config["test_predictions"] = str(ROOT / "predictions/test_predictions.csv")
config["report"] = str(report_path)
config_path.write_text(json.dumps(config, indent=2, allow_nan=False), encoding="utf-8")
print(report_path)
# END REGISTERED SOURCE BLOCK


#### Earlier methodology setup (cell 1)

In [104]:
%%project_source historical/v2/methodology_gap_analysis_v2.ipynb::cell1 0
from pathlib import Path
import json, hashlib, math, warnings
import numpy as np
import pandas as pd
import matplotlib.pyplot as plt
from PIL import Image
from scipy.fft import dctn
from scipy.stats import chi2_contingency
from sklearn.calibration import calibration_curve
from sklearn.linear_model import LogisticRegression
from sklearn.metrics import (
    accuracy_score, precision_score, recall_score, f1_score,
    roc_auc_score, average_precision_score, brier_score_loss,
    log_loss, confusion_matrix
)
from sklearn.model_selection import train_test_split

ORIGINAL_ROOT = Path(r"F:\data sci\project\multimodal-fake-news-detection").resolve()
V2_ROOT = Path(r"F:\data sci\project\v2").resolve()
OUTPUT_ROOT = V2_ROOT / "outputs"
MANIFEST_ROOT = V2_ROOT / "manifests"
RAW_ROOT = ORIGINAL_ROOT / "data" / "raw" / "fakeddit"
PROCESSED_ROOT = ORIGINAL_ROOT / "data" / "processed" / "fakeddit"
RESULTS_ROOT = ORIGINAL_ROOT / "results"
SEED = 2026

assert ORIGINAL_ROOT.exists(), ORIGINAL_ROOT
assert V2_ROOT != ORIGINAL_ROOT and ORIGINAL_ROOT not in V2_ROOT.parents
OUTPUT_ROOT.mkdir(parents=True, exist_ok=True)
MANIFEST_ROOT.mkdir(parents=True, exist_ok=True)

def save_json(name, obj):
    path = OUTPUT_ROOT / name
    path.write_text(json.dumps(obj, indent=2, default=str), encoding="utf-8")
    return path

def raw_path(split):
    name = {"train":"multimodal_train.tsv", "validation":"multimodal_validate.tsv", "test":"multimodal_test_public.tsv"}[split]
    return RAW_ROOT / "multimodal_only_samples" / name

def read_raw(split, columns=None):
    return pd.read_csv(raw_path(split), sep="\t", usecols=columns, low_memory=False)

def metrics(y, p, threshold=0.5):
    y = np.asarray(y, dtype=int); p = np.clip(np.asarray(p, dtype=float), 1e-7, 1-1e-7)
    pred = (p >= threshold).astype(int)
    return {
        "n": int(len(y)), "threshold": float(threshold),
        "accuracy": float(accuracy_score(y, pred)),
        "precision": float(precision_score(y, pred, zero_division=0)),
        "recall": float(recall_score(y, pred, zero_division=0)),
        "f1": float(f1_score(y, pred, zero_division=0)),
        "macro_f1": float(f1_score(y, pred, average="macro", zero_division=0)),
        "roc_auc": float(roc_auc_score(y, p)) if len(np.unique(y)) == 2 else np.nan,
        "pr_auc": float(average_precision_score(y, p)) if len(np.unique(y)) == 2 else np.nan,
        "brier": float(brier_score_loss(y, p)),
        "log_loss": float(log_loss(y, p, labels=[0,1])),
        "confusion_matrix": confusion_matrix(y, pred, labels=[0,1]).tolist(),
    }

print("Original (read-only):", ORIGINAL_ROOT)
print("v2 outputs:", V2_ROOT)
# END REGISTERED SOURCE BLOCK


### Recorded configuration and dependencies

These are recorded project settings and environment snapshots, not a promise that every pinned version installs on every platform. Use a compatible Python/PyTorch/torchvision environment for the available hardware. The ordinary and source-disjoint configurations belong to different experiments.

#### `multimodal-fake-news-detection/configs/base.yaml`

```
project:
  name: multimodal-fake-news-detection
  seed: 42

task:
  type: binary_classification
  num_classes: 2

data:
  train_ratio: 0.70
  validation_ratio: 0.15
  test_ratio: 0.15
  num_workers: 4

training:
  epochs: 5
  early_stopping_patience: 2

evaluation:
  metrics:
    - accuracy
    - precision
    - recall
    - f1
    - roc_auc
    - pr_auc

```

#### `multimodal-fake-news-detection/configs/fakeddit_data.yaml`

```
dataset:
  name: fakeddit
  version: "2.0"
  task: binary_classification
  source_label_column: 2_way_label

development_subset:
  seed: 42

  original:
    train: 20000
    validation: 3000
    test: 3000

  cleaned_multimodal:
    train: 13129
    validation: 1962
    test: 1965

paths:
  train: data/processed/fakeddit/development_clean/train.parquet
  validation: data/processed/fakeddit/development_clean/validation.parquet
  test: data/processed/fakeddit/development_clean/test.parquet

modalities:
  text:
    column: text
    source: clean_title

  image:
    column: image_path
    root: data/raw/fakeddit/development_images

cleaning:
  require_existing_image: true
  require_valid_image: true

  excluded_placeholder:
    sha256: faa24ec881e6040655c187a681d6dc496eb8aa41e1bd0652a180b3a40b457187
    source_subreddit: psbattle_artwork
    reason: repeated regional-unavailable placeholder image

splits:
  preserve_official_fakeddit_boundaries: true
  identical_sample_ids_across_modalities: true

text_processing:
  tokenizer: roberta-base
  max_length: 64

evaluation:
  main_metrics:
    - accuracy
    - precision
    - recall
    - f1
    - roc_auc
    - pr_auc

notes:
  class_distribution_shift_after_image_filtering: true
  placeholder_images_are_class_conditional: true
  do_not_rebalance_main_benchmark: true

```

#### `multimodal-fake-news-detection/requirements.txt`

```
accelerate==1.14.0
aiohappyeyeballs==2.7.1
aiohttp==3.14.3
aiosignal==1.4.0
annotated-doc==0.0.5
anyio==4.14.2
argon2-cffi==25.1.0
argon2-cffi-bindings==26.1.0
arrow==1.4.0
asttokens==3.0.2
async-lru==2.3.0
attrs==26.1.0
babel==2.18.0
beautifulsoup4==4.15.0
bleach==6.4.0
certifi==2026.7.22
cffi==2.1.1
charset-normalizer==3.5.1
click==8.5.0
cloudpickle==3.1.2
colorama==0.4.6
comm==0.2.3
contourpy==1.3.3
cycler==0.12.1
datasets==5.0.1
debugpy==1.8.21
defusedxml==0.7.1
dill==0.4.1
executing==2.2.1
fastjsonschema==2.22.2
filelock==3.32.5
fonttools==4.64.0
fqdn==1.5.1
frozenlist==1.8.0
fsspec==2026.6.0
gdown==6.1.0
h11==0.16.0
hf-xet==1.6.0
httpcore==1.0.9
httpx==0.28.1
huggingface_hub==1.29.0
idna==3.19
iniconfig==2.3.0
ipykernel==7.3.0
ipython==9.17.0
ipython_pygments_lexers==1.1.1
isoduration==20.11.0
jedi==0.20.0
Jinja2==3.1.6
joblib==1.6.0
json5==0.15.0
jsonpointer==3.1.1
jsonschema==4.26.0
jsonschema-specifications==2025.9.1
jupyter-events==0.12.1
jupyter-lsp==2.3.1
jupyter_builder==1.2.2
jupyter_client==8.10.0
jupyter_core==5.9.1
jupyter_server==2.21.0
jupyter_server_terminals==0.5.4
jupyterlab==4.6.3
jupyterlab_pygments==0.3.0
jupyterlab_server==2.28.0
kiwisolver==1.5.1
lark==1.3.1
lightning-utilities==0.15.3
markdown-it-py==4.2.0
MarkupSafe==3.0.3
matplotlib==3.11.1
matplotlib-inline==0.2.2
mdurl==0.1.2
mistune==3.3.4
mpmath==1.3.0
multidict==6.7.1
multiprocess==0.70.19
narwhals==2.25.0
nbclient==0.11.0
nbconvert==7.17.1
nbformat==5.11.1
nest-asyncio2==1.7.2
networkx==3.6.1
notebook_shim==0.2.4
numpy==2.5.2
opencv-python==5.0.0.93
packaging==26.3
pandas==3.0.5
pandocfilters==1.5.1
parso==0.8.7
pillow==12.3.0
platformdirs==4.11.5
pluggy==1.6.0
prometheus_client==0.26.0
prompt_toolkit==3.0.53
propcache==0.5.2
psutil==7.2.2
pure_eval==0.2.3
pyarrow==25.0.1
pycparser==3.0
Pygments==2.21.0
pyparsing==3.3.2
PySocks==1.7.1
pytest==9.1.1
python-dateutil==2.9.0.post0
python-dotenv==1.2.3
python-json-logger==4.2.0
pywinpty==3.0.5
PyYAML==6.0.3
pyzmq==27.2.0
referencing==0.37.0
regex==2026.8.31
requests==2.34.2
rfc3339-validator==0.1.4
rfc3986-validator==0.1.1
rfc3987-syntax==1.1.0
rich==15.0.0
rpds-py==2026.6.3
safetensors==0.8.0
scikit-learn==1.9.0
scipy==1.18.1
Send2Trash==2.1.0
setuptools==84.0.0
shellingham==1.5.4
six==1.17.0
soupsieve==2.9.2
stack-data==0.6.3
sympy==1.14.0
terminado==0.18.1
threadpoolctl==3.6.0
timm==1.0.29
tinycss2==1.5.1
tokenizers==0.23.1
torch==2.13.0
torchaudio==2.11.0
torchmetrics==1.9.0
torchvision==0.28.0
tornado==6.5.8
tqdm==4.70.0
traitlets==5.16.1
transformers==5.16.1
typer==0.27.2
typing_extensions==4.16.0
tzdata==2026.3
uri-template==1.3.0
urllib3==2.7.0
wcwidth==0.8.3
webcolors==25.10.0
webencodings==0.6.1
websocket-client==1.9.2
xxhash==4.0.1
yarl==1.24.5

```

#### `multimodal-fake-news-detection/requirements-desktop.txt`

```
accelerate==1.14.0
aiohappyeyeballs==2.7.1
aiohttp==3.14.3
aiosignal==1.4.0
annotated-doc==0.0.5
anyio==4.14.2
argon2-cffi==25.1.0
argon2-cffi-bindings==26.1.0
arrow==1.4.0
asttokens==3.0.2
async-lru==2.3.0
attrs==26.1.0
babel==2.18.0
beautifulsoup4==4.15.0
bleach==6.4.0
certifi==2026.7.22
cffi==2.1.1
charset-normalizer==3.5.1
click==8.5.0
cloudpickle==3.1.2
colorama==0.4.6
comm==0.2.3
contourpy==1.3.3
cycler==0.12.1
datasets==5.0.1
debugpy==1.8.21
defusedxml==0.7.1
dill==0.4.1
executing==2.2.1
fastjsonschema==2.22.2
filelock==3.32.5
fonttools==4.64.0
fqdn==1.5.1
frozenlist==1.8.0
fsspec==2026.6.0
gdown==6.1.0
h11==0.16.0
hf-xet==1.6.0
httpcore==1.0.9
httpx==0.28.1
huggingface_hub==1.29.0
idna==3.19
iniconfig==2.3.0
ipykernel==7.3.0
ipython==9.17.0
ipython_pygments_lexers==1.1.1
isoduration==20.11.0
jedi==0.20.0
Jinja2==3.1.6
joblib==1.6.0
json5==0.15.0
jsonpointer==3.1.1
jsonschema==4.26.0
jsonschema-specifications==2025.9.1
jupyter-events==0.12.1
jupyter-lsp==2.3.1
jupyter_builder==1.2.2
jupyter_client==8.10.0
jupyter_core==5.9.1
jupyter_server==2.21.0
jupyter_server_terminals==0.5.4
jupyterlab==4.6.3
jupyterlab_pygments==0.3.0
jupyterlab_server==2.28.0
kiwisolver==1.5.1
lark==1.3.1
lightning-utilities==0.15.3
markdown-it-py==4.2.0
MarkupSafe==3.0.3
matplotlib==3.11.1
matplotlib-inline==0.2.2
mdurl==0.1.2
mistune==3.3.4
mpmath==1.3.0
multidict==6.7.1
multiprocess==0.70.19
narwhals==2.25.0
nbclient==0.11.0
nbconvert==7.17.1
nbformat==5.11.1
nest-asyncio2==1.7.2
networkx==3.6.1
notebook_shim==0.2.4
numpy==2.5.2
opencv-python==5.0.0.93
packaging==26.3
pandas==3.0.5
pandocfilters==1.5.1
parso==0.8.7
pillow==12.3.0
platformdirs==4.11.5
pluggy==1.6.0
prometheus_client==0.26.0
prompt_toolkit==3.0.53
propcache==0.5.2
psutil==7.2.2
pure_eval==0.2.3
pyarrow==25.0.1
pycparser==3.0
Pygments==2.21.0
pyparsing==3.3.2
PySocks==1.7.1
pytest==9.1.1
python-dateutil==2.9.0.post0
python-dotenv==1.2.3
python-json-logger==4.2.0
pywinpty==3.0.5
PyYAML==6.0.3
pyzmq==27.2.0
referencing==0.37.0
regex==2026.8.31
requests==2.34.2
rfc3339-validator==0.1.4
rfc3986-validator==0.1.1
rfc3987-syntax==1.1.0
rich==15.0.0
rpds-py==2026.6.3
safetensors==0.8.0
scikit-learn==1.9.0
scipy==1.18.1
Send2Trash==2.1.0
setuptools==84.0.0
shellingham==1.5.4
six==1.17.0
soupsieve==2.9.2
stack-data==0.6.3
sympy==1.14.0
terminado==0.18.1
threadpoolctl==3.6.0
timm==1.0.29
tinycss2==1.5.1
tokenizers==0.23.1
torchmetrics==1.9.0
tornado==6.5.8
tqdm==4.70.0
traitlets==5.16.1
transformers==5.16.1
typer==0.27.2
typing_extensions==4.16.0
tzdata==2026.3
uri-template==1.3.0
urllib3==2.7.0
wcwidth==0.8.3
webcolors==25.10.0
webencodings==0.6.1
websocket-client==1.9.2
xxhash==4.0.1
yarl==1.24.5

```

#### `v2/experiments/source_disjoint/experiment_config.json`

```
{
  "experiment": "source_disjoint",
  "created_utc": "2026-09-15T11:18:00.664633+00:00",
  "seed": 42,
  "project_root": "F:\\data sci\\project\\multimodal-fake-news-detection",
  "source_manifest": "F:\\data sci\\project\\v2\\manifests\\source_disjoint.parquet",
  "isolated_manifest": "F:\\data sci\\project\\v2\\experiments\\source_disjoint\\manifests\\source_disjoint.parquet",
  "manifest_sha256": "f7feb3531ef6decd1ea95af9dce8eeb7dbf7d2f7670b8db68c614a721308cc52",
  "split_counts": {
    "train": 10524,
    "validation": 3793,
    "test": 2739
  },
  "positive_class": 1,
  "classification_threshold": 0.5,
  "roberta": {
    "base_model": "roberta-base",
    "pretrained_base_weights": true,
    "max_length": 64,
    "batch_size": 16,
    "optimizer": "AdamW",
    "learning_rate": 2e-05,
    "weight_decay": 0.01,
    "gradient_clipping": 1.0,
    "warmup_fraction": 0.1,
    "max_epochs": 3,
    "selection_metric": "validation_macro_f1",
    "checkpoint": "F:\\data sci\\project\\v2\\experiments\\source_disjoint\\checkpoints\\roberta"
  },
  "resnet50": {
    "base_model": "resnet50",
    "weights": "IMAGENET1K_V2",
    "fine_tune": "full network",
    "input_size": [
      224,
      224
    ],
    "batch_size": 32,
    "optimizer": "AdamW",
    "learning_rate": 0.0001,
    "weight_decay": 0.01,
    "max_epochs": 3,
    "selection_metric": "validation_macro_f1",
    "checkpoint": "F:\\data sci\\project\\v2\\experiments\\source_disjoint\\checkpoints\\resnet50\\best_model.pt"
  },
  "fusion": {
    "formula": "alpha * p_text + (1 - alpha) * p_image",
    "alpha_search": [
      0.0,
      0.05,
      0.1,
      0.15,
      0.2,
      0.25,
      0.3,
      0.35,
      0.4,
      0.45,
      0.5,
      0.55,
      0.6,
      0.65,
      0.7,
      0.75,
      0.8,
      0.85,
      0.9,
      0.95,
      1.0
    ],
    "selection_metric": "validation_macro_f1",
    "tie_break": "closest to 0.50, then lower alpha",
    "selected_alpha": 0.0,
    "locked_utc": "2026-09-15T11:28:39.694083+00:00"
  },
  "calibration": {
    "ece_bins": 10,
    "convention": "confidence bins from 0.5 to 1.0"
  },
  "bootstrap": {
    "iterations": 5000,
    "seed": 42,
    "paired": true
  },
  "packages": {
    "python": "3.12.3",
    "torch": "2.13.0+cu126",
    "torchvision": "0.28.0+cu126",
    "transformers": "5.16.1",
    "pandas": "3.0.5",
    "numpy": "2.5.2",
    "scikit_learn": "1.9.0",
    "scipy": "1.18.1"
  },
  "hardware": {
    "cuda_available": true,
    "cuda_version": "12.6",
    "gpu": "NVIDIA GeForce RTX 2070 SUPER"
  },
  "test_evaluated_utc": "2026-09-15T11:33:30.919858+00:00",
  "test_predictions": "F:\\data sci\\project\\v2\\experiments\\source_disjoint\\predictions\\test_predictions.csv",
  "report": "F:\\data sci\\project\\v2\\experiments\\source_disjoint\\reports\\source_disjoint_results.md"
}
```

<a id="reproduce"></a>
## 11. Saved evidence and reproduction controls

The next collapsed cell stores a compressed copy of the saved evidence, including predictions and manifests. It is data, not a trained model or hidden implementation. All Python implementation is visible above. The archive is extracted only into a fresh directory, and filenames are checked before extraction. No original project file is modified.

In [105]:
EVIDENCE_ARCHIVE_B64 = '...'
EXPECTED_SOURCE_HASHES = {'multimodal-fake-news-detection/scripts/audit_fakeddit.py': 'd4fd48d8cc076a2452dd35607d77bf6a57ead41491d7f6371ea57186b0d551a7', 'multimodal-fake-news-detection/scripts/audit_split_leakage.py': '47fe810833df421065be9ea249c68b5741608780fefd7c5fb90b2e0f75ff52b9', 'multimodal-fake-news-detection/scripts/prepare_fakeddit.py': 'be2a99e0a7ba9378453bbeebe4db45e2f80573fc58cec88fc2927e81b1b634c4', 'multimodal-fake-news-detection/scripts/create_dev_subset.py': '83d207a45502c8fa5196fa80bd0a645833cec1b0f61051ecec914c55cb4a3557', 'multimodal-fake-news-detection/scripts/download_dev_images.py': '03b09707f152859b110a5772994866d744adc3a43e1a19137727e7ef5941fa57', 'multimodal-fake-news-detection/scripts/audit_image_integrity.py': '023e7d1d1db932c160fb5718df72e893209c4a0495a74ba89d5e99d6776cd0cf', 'multimodal-fake-news-detection/scripts/inspect_duplicate_hashes.py': 'bf92a068c85a216817f098ba9ae072012117d822899700fe06be587b97373ca7', 'multimodal-fake-news-detection/scripts/create_clean_multimodal_manifests.py': 'f197933f57c4c730b0fab509c145d655afd1c018f854b23e07a22b969111645a', 'multimodal-fake-news-detection/scripts/analyse_placeholder_sources.py': '2a3ea9df3e7e85bb6bbf6ad21e9c5545ea2f1c1aa374eb0560f3154f9e33a57f', 'multimodal-fake-news-detection/scripts/freeze_fakeddit_data.py': 'e28103c32e39fdc972d2e767503455b5ce438ea70da0e1463b156b0c612ea154', 'multimodal-fake-news-detection/scripts/generate_eda_figures.py': '3f70f7b5dfa8ee16ab892c3f900f8f4d69e6536dcb0cf19dd3e10beaad0071a5', 'multimodal-fake-news-detection/scripts/audit_token_lengths.py': '6804b08ffafea755f52c6c126e7a5dab0495b86d927221dfd60e10ce75526799', 'multimodal-fake-news-detection/scripts/train_roberta_baseline.py': '13684f20c54175060ea306d60641f065000dc1ce61ae18e1a0e95e1973906091', 'multimodal-fake-news-detection/scripts/plot_roberta_baseline.py': '96d9e87cc106fdefcdf9b2548c7c86c8153d333e5940aea9e288c3d02cfef202', 'multimodal-fake-news-detection/scripts/train_resnet_baseline.py': 'a8f7e21493c7d391b6c3013ee1212054b1bd590cf5fc8b47a9ce99293d988f8f', 'multimodal-fake-news-detection/scripts/extract_multimodal_features.py': 'f9fbcc5f6ccbedcb7e8c7064bcfd17de48a89582537851dafdbc3e54504cb665', 'multimodal-fake-news-detection/scripts/train_multimodal_fusion.py': '3e68497230c7e422e4cad06e513b4ea38843554d01e99a4ea9cf47b7e6f881e3', 'multimodal-fake-news-detection/scripts/tune_multimodal_fusion.py': 'd43899356ca268691114683c6c7dd7a2d0d2903915005d9457c70a110d3ff7bd', 'multimodal-fake-news-detection/scripts/evaluate_linear_fusion.py': '0738418c3c8befe5a8fb932a3eb220be58d8d8390f84d29f5967f17928da6ec7', 'multimodal-fake-news-detection/scripts/export_baseline_probabilities.py': 'a89f4a953b215ad1a30a38bd612f29fde83ec24ef3789fcbd4e2f3cd3f52bf99', 'multimodal-fake-news-detection/scripts/evaluate_late_fusion.py': 'afd48c5d789e045a1d918e89e0f91061cf71197a341efbb56a792d39a5f9017f', 'multimodal-fake-news-detection/scripts/compare_fusion_vs_roberta.py': '9d45a57e1a997c14ce4e5ee8dd5394b52835e07ac7a4dec42db886103e68a07f', 'multimodal-fake-news-detection/scripts/analyse_calibration.py': '7f2a89322f5adfad2d0687751673d710c54eca1632e2c5da38223eba4b1556ed', 'multimodal-fake-news-detection/scripts/analyse_missing_modality.py': '2f733b24d2560a5b398e6b50b1d6f7254192d93c02837ab7b0fb724b17ec9dd7', 'multimodal-fake-news-detection/scripts/analyse_model_errors.py': '9b07320810e0f0ac93f8d49b4a6414902f70781501d09fd515605410d42e7988', 'multimodal-fake-news-detection/scripts/generate_roberta_shap_cases.py': '175303ca5e803ad1575fdf628226006fb0d164ace87206877347bfca21e1a171', 'multimodal-fake-news-detection/scripts/generate_gradcam_cases.py': 'e3b2285679cb0e1063d5916362ecd290382017b2699a9f4f9b9a77d6439b0524', 'multimodal-fake-news-detection/scripts/build_multimodal_case_studies.py': '80798863bd55b16a1b2619bf0486ef118e66936d9f7c7f954f46511b30d17933', 'multimodal-fake-news-detection/scripts/create_final_holdout_candidates.py': '6680ea2826211949f1eb28e1e7ebc0d8c0748abc2986e36e7ea5cd4a8c039cec', 'multimodal-fake-news-detection/scripts/prepare_final_holdout.py': '7d358b12eb6d4a657a75818f62469347d0b1f0d80a1b14ea6ae7d2572fbd05d6', 'multimodal-fake-news-detection/scripts/evaluate_final_holdout.py': 'f840fad628de5b07152e4dec74790045dacdd1881d03e2e96d8b62112f33b83f', 'v2/methodology_gap_analysis_v2.ipynb::cell1': 'd0e55062350d96b01db14aeef14edf258760be54b28a64b9d530037d0331f40f', 'v2/methodology_gap_analysis_v2.ipynb::cell3': '47f157225242fe0c83da57eb9b9f671501ff675e686845ac82bbdea96a6c0be3', 'v2/methodology_gap_analysis_v2.ipynb::cell5': 'a311a9a7725d11b02bcf7d66630efc49881f487f09269691dbaf89cdbad6ec6d', 'v2/methodology_gap_analysis_v2.ipynb::cell7': 'e3c611fe46fa0558a751959e1a3ca5016315d25d91727abee5214ad17fd2d988', 'v2/methodology_gap_analysis_v2.ipynb::cell9': '5d0d21664e7a44cdb0356c3b04220e6aa1417f911edd7721c106cf29e5023db6', 'v2/methodology_gap_analysis_v2.ipynb::cell11': '7ea08042e1e81898d9325b6077be12983da73961f4a1c2b2f2f4682992b052aa', 'v2/methodology_gap_analysis_v2.ipynb::cell13': '636fe14733ece2e26ccb781d38c014ac803b9c5ee06c2752d7ad5e2110ef2bc6', 'v2/methodology_gap_analysis_v2.ipynb::cell15': 'df75c7bf8f664768f06713353924656b7b5e2e164aac0c829888b1faea176c53', 'v2/experiments/source_disjoint/run_source_disjoint.py': 'daa0441868b2c7c565ac0053813809c2dcd1e708ca2d7a4a6097a82f00f57388', 'tools/verify_saved_results.py': 'ce1b28e97eadba802c58130084962d78eaa4f9262f8f240773b533dff2a6cf6e', 'multimodal-fake-news-detection/tests/test_environment.py': '58e03bfdda67d360be291ffebc885383ee597da22d2e856ceb93a96031d1a033', 'multimodal-fake-news-detection/src/fake_news/__init__.py': '01ba4719c80b6fe911b091a7c05124b64eeece964e09c058ef8f9805daca546b', 'multimodal-fake-news-detection/src/fake_news/data/__init__.py': '01ba4719c80b6fe911b091a7c05124b64eeece964e09c058ef8f9805daca546b', 'multimodal-fake-news-detection/src/fake_news/evaluation/__init__.py': '01ba4719c80b6fe911b091a7c05124b64eeece964e09c058ef8f9805daca546b', 'multimodal-fake-news-detection/src/fake_news/explainability/__init__.py': '01ba4719c80b6fe911b091a7c05124b64eeece964e09c058ef8f9805daca546b', 'multimodal-fake-news-detection/src/fake_news/models/__init__.py': '01ba4719c80b6fe911b091a7c05124b64eeece964e09c058ef8f9805daca546b', 'multimodal-fake-news-detection/src/fake_news/training/__init__.py': '01ba4719c80b6fe911b091a7c05124b64eeece964e09c058ef8f9805daca546b', 'historical/v2/experiments/source_disjoint/run_source_disjoint.py': '36acc2b421bd831702cb09d4293e12f6090c21e522a3290b82031fb253c7caad', 'historical/v2/experiments/source_disjoint/build_report.py': '11d3641acc8886bdadfaa2d24e480b4ebfac5388f7140e112d6f07107a534468', 'historical/v2/methodology_gap_analysis_v2.ipynb::cell1': 'b20975653e1232fc2e592046405f541f00b11b8a4025723996388811038087fd'}
NOTEBOOK_DOCUMENTS = {'v2/methodology_gap_analysis_v2.ipynb': {'cells': [{'cell_type': 'markdown', 'id': '4e390fca', 'metadata': {}, 'source': ['# Fakeddit multimodal methodology audit — v2\n', '\n', 'This notebook adds the methodological checks that were missing from the original project while preserving the original code, data, checkpoints, and results. It reads from the sibling `multimodal-fake-news-detection` folder and writes only to this `v2` folder.\n', '\n', 'The notebook covers:\n', '\n', '1. binary-label semantics and internal consistency;\n', '2. class-dependent image-selection bias;\n', '3. a fairer validation-tuned and calibrated RoBERTa comparison;\n', '4. source, domain, and time subgroup performance plus a source-only shortcut baseline;\n', '5. perceptual-image duplicate screening;\n', '6. source-disjoint and chronological manifests for stronger future retraining;\n', '7. explainability coverage and reporting consistency checks.\n', '\n', 'The final holdout is used only for locked evaluation of predeclared controls. No original model or result is overwritten.']}, {'cell_type': 'code', 'execution_count': None, 'id': '150aecf6', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:48.042916Z', 'iopub.status.busy': '2026-09-09T12:46:48.041916Z', 'iopub.status.idle': '2026-09-09T12:46:49.845246Z', 'shell.execute_reply': '2026-09-09T12:46:49.845246Z'}}, 'outputs': [], 'source': ['from pathlib import Path\n', 'import json, hashlib, math, warnings\n', 'import numpy as np\n', 'import pandas as pd\n', 'import matplotlib.pyplot as plt\n', 'from PIL import Image\n', 'from scipy.fft import dctn\n', 'from scipy.stats import chi2_contingency\n', 'from sklearn.calibration import calibration_curve\n', 'from sklearn.linear_model import LogisticRegression\n', 'from sklearn.metrics import (\n', '    accuracy_score, precision_score, recall_score, f1_score,\n', '    roc_auc_score, average_precision_score, brier_score_loss,\n', '    log_loss, confusion_matrix\n', ')\n', 'from sklearn.model_selection import train_test_split\n', '\n', '# Open the notebook from v2 or the submission repository root.\n', 'REPO_ROOT = Path.cwd().resolve()\n', 'if REPO_ROOT.name == "v2":\n', '    REPO_ROOT = REPO_ROOT.parent\n', 'ORIGINAL_ROOT = REPO_ROOT / "multimodal-fake-news-detection"\n', 'V2_ROOT = REPO_ROOT / "v2"\n', 'OUTPUT_ROOT = V2_ROOT / "outputs"\n', 'MANIFEST_ROOT = V2_ROOT / "manifests"\n', 'RAW_ROOT = ORIGINAL_ROOT / "data" / "raw" / "fakeddit"\n', 'PROCESSED_ROOT = ORIGINAL_ROOT / "data" / "processed" / "fakeddit"\n', 'RESULTS_ROOT = ORIGINAL_ROOT / "results"\n', 'SEED = 2026\n', '\n', 'assert ORIGINAL_ROOT.exists(), ORIGINAL_ROOT\n', 'assert V2_ROOT != ORIGINAL_ROOT and ORIGINAL_ROOT not in V2_ROOT.parents\n', 'OUTPUT_ROOT.mkdir(parents=True, exist_ok=True)\n', 'MANIFEST_ROOT.mkdir(parents=True, exist_ok=True)\n', '\n', 'def save_json(name, obj):\n', '    path = OUTPUT_ROOT / name\n', '    path.write_text(json.dumps(obj, indent=2, default=str), encoding="utf-8")\n', '    return path\n', '\n', 'def raw_path(split):\n', '    name = {"train":"multimodal_train.tsv", "validation":"multimodal_validate.tsv", "test":"multimodal_test_public.tsv"}[split]\n', '    return RAW_ROOT / "multimodal_only_samples" / name\n', '\n', 'def read_raw(split, columns=None):\n', '    return pd.read_csv(raw_path(split), sep="\\t", usecols=columns, low_memory=False)\n', '\n', 'def metrics(y, p, threshold=0.5):\n', '    y = np.asarray(y, dtype=int); p = np.clip(np.asarray(p, dtype=float), 1e-7, 1-1e-7)\n', '    pred = (p >= threshold).astype(int)\n', '    return {\n', '        "n": int(len(y)), "threshold": float(threshold),\n', '        "accuracy": float(accuracy_score(y, pred)),\n', '        "precision": float(precision_score(y, pred, zero_division=0)),\n', '        "recall": float(recall_score(y, pred, zero_division=0)),\n', '        "f1": float(f1_score(y, pred, zero_division=0)),\n', '        "macro_f1": float(f1_score(y, pred, average="macro", zero_division=0)),\n', '        "roc_auc": float(roc_auc_score(y, p)) if len(np.unique(y)) == 2 else np.nan,\n', '        "pr_auc": float(average_precision_score(y, p)) if len(np.unique(y)) == 2 else np.nan,\n', '        "brier": float(brier_score_loss(y, p)),\n', '        "log_loss": float(log_loss(y, p, labels=[0,1])),\n', '        "confusion_matrix": confusion_matrix(y, pred, labels=[0,1]).tolist(),\n', '    }\n', '\n', 'print("Original (read-only):", ORIGINAL_ROOT)\n', 'print("v2 outputs:", V2_ROOT)']}, {'cell_type': 'markdown', 'id': '4d875460', 'metadata': {}, 'source': ['## 1. Verify label semantics\n', '\n', "Fakeddit's six-way label `0` is the true-content category; the other five categories are forms of false or misleading content. The binary encoding is therefore checked programmatically: binary class `1` must correspond exactly to six-way class `0`, and binary class `0` to six-way classes `1–5`."]}, {'cell_type': 'code', 'execution_count': None, 'id': 'cf69b2b5', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:49.847787Z', 'iopub.status.busy': '2026-09-09T12:46:49.846782Z', 'iopub.status.idle': '2026-09-09T12:46:51.906215Z', 'shell.execute_reply': '2026-09-09T12:46:51.906215Z'}}, 'outputs': [], 'source': ['label_rows = []\n', 'label_tables = {}\n', 'for split in ["train", "validation", "test"]:\n', '    d = read_raw(split, ["id", "2_way_label", "3_way_label", "6_way_label"])\n', '    tab = pd.crosstab(d["2_way_label"], d["6_way_label"])\n', '    label_tables[split] = tab\n', '    consistent = ((d["2_way_label"] == 1) == (d["6_way_label"] == 0))\n', '    label_rows.append({\n', '        "split": split, "n": len(d), "consistent_n": int(consistent.sum()),\n', '        "inconsistent_n": int((~consistent).sum()), "consistent_pct": float(100*consistent.mean())\n', '    })\n', '    display(tab)\n', '\n', 'label_audit = pd.DataFrame(label_rows)\n', 'label_audit.to_csv(OUTPUT_ROOT / "label_semantics_audit.csv", index=False)\n', 'assert label_audit["inconsistent_n"].sum() == 0\n', 'semantics = {\n', '    "binary_class_1": "true/real content",\n', '    "binary_class_0": "fake or misleading content (six-way classes 1-5)",\n', '    "verification": label_rows,\n', '    "limitation": "This verifies dataset encoding, not the factual correctness of every distant-supervision label."\n', '}\n', 'save_json("label_semantics.json", semantics)\n', 'display(label_audit)']}, {'cell_type': 'markdown', 'id': '3a8ba1ee', 'metadata': {}, 'source': ['## 2. Quantify selection bias caused by image availability\n', '\n', 'Equal sample IDs make comparisons between modalities fair within the retained subset. They do not make that subset representative. This section measures retention by label, year, domain, and subreddit and tests whether retention is independent of the binary label.']}, {'cell_type': 'code', 'execution_count': None, 'id': 'de8fac17', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:51.908257Z', 'iopub.status.busy': '2026-09-09T12:46:51.908257Z', 'iopub.status.idle': '2026-09-09T12:46:55.460716Z', 'shell.execute_reply': '2026-09-09T12:46:55.460716Z'}}, 'outputs': [], 'source': ['status_parts = []\n', 'for split in ["train", "validation", "test"]:\n', '    p = PROCESSED_ROOT / "development_clean" / f"{split}_with_image_status.parquet"\n', '    s = pd.read_parquet(p)\n', '    meta = read_raw(split, ["id", "subreddit", "domain", "created_utc", "2_way_label"])\n', '    s["id"] = s["id"].astype(str); meta["id"] = meta["id"].astype(str)\n', '    s = s.merge(meta, on="id", how="left", validate="one_to_one")\n', '    s["retained"] = s["image_usable"].fillna(False).astype(bool)\n', '    s["year"] = pd.to_datetime(s["created_utc"], unit="s", errors="coerce", utc=True).dt.year\n', '    status_parts.append(s)\n', 'status = pd.concat(status_parts, ignore_index=True)\n', '\n', 'retention = (status.groupby(["split", "label"])["retained"]\n', '             .agg(total="size", retained="sum", retention_rate="mean").reset_index())\n', 'retention["removed"] = retention["total"] - retention["retained"]\n', 'retention.to_csv(OUTPUT_ROOT / "selection_retention_by_label.csv", index=False)\n', '\n', 'contingency = pd.crosstab(status["label"], status["retained"])\n', 'chi2, p_value, _, _ = chi2_contingency(contingency)\n', 'n = contingency.to_numpy().sum()\n', 'cramers_v = math.sqrt(chi2 / n)\n', 'bias_summary = {\n', '    "n": int(n), "chi_square": float(chi2), "p_value": float(p_value),\n', '    "cramers_v": float(cramers_v),\n', '    "interpretation": "Large dependence means complete-case filtering changes the target population. Macro-F1 does not remove this selection bias."\n', '}\n', 'save_json("selection_bias_summary.json", bias_summary)\n', '\n', 'for group in ["subreddit", "domain", "year"]:\n', '    g = (status.groupby(group, dropna=False)["retained"]\n', '         .agg(total="size", retained="sum", retention_rate="mean").reset_index())\n', '    g["removed"] = g["total"] - g["retained"]\n', '    g.sort_values(["total", "retention_rate"], ascending=[False, True]).to_csv(\n', '        OUTPUT_ROOT / f"selection_retention_by_{group}.csv", index=False)\n', '\n', 'display(retention)\n', 'print(bias_summary)\n', '\n', 'fig, ax = plt.subplots(figsize=(7,4))\n', 'for split, grp in retention.groupby("split"):\n', '    ax.plot(grp["label"].astype(str), grp["retention_rate"], marker="o", label=split)\n', 'ax.set(xlabel="Binary label (0=fake/misleading, 1=true)", ylabel="Image retention rate", ylim=(0,1),\n', '       title="Image filtering is strongly class-dependent")\n', 'ax.legend(); fig.tight_layout()\n', 'fig.savefig(OUTPUT_ROOT / "selection_retention_by_label.png", dpi=180)\n', 'plt.show()']}, {'cell_type': 'markdown', 'id': '0e54206c', 'metadata': {}, 'source': ['## 3. Fair text-only threshold and calibration controls\n', '\n', 'The original fusion weight was selected on validation macro-F1 while RoBERTa used the default 0.5 threshold. This section gives RoBERTa the same opportunity to tune its decision threshold. It also fits Platt calibration on one stratified half of validation and selects its threshold on the other half, then evaluates each predeclared variant once on the frozen holdout.']}, {'cell_type': 'code', 'execution_count': None, 'id': '6fe2166a', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:55.462761Z', 'iopub.status.busy': '2026-09-09T12:46:55.462761Z', 'iopub.status.idle': '2026-09-09T12:46:58.608870Z', 'shell.execute_reply': '2026-09-09T12:46:58.608870Z'}}, 'outputs': [], 'source': ['val = pd.read_csv(RESULTS_ROOT / "metrics" / "baseline_probabilities" / "roberta_validation.csv")\n', 'final = pd.read_csv(RESULTS_ROOT / "metrics" / "final_evaluation" / "final_predictions.csv")\n', 'val = val.rename(columns={"probability_class_1":"p_text"})\n', '\n', 'threshold_grid = np.linspace(0.05, 0.95, 181)\n', 'threshold_scores = pd.DataFrame({\n', '    "threshold": threshold_grid,\n', '    "validation_macro_f1": [metrics(val.label, val.p_text, t)["macro_f1"] for t in threshold_grid]\n', '})\n', 'best_t = float(threshold_scores.sort_values(["validation_macro_f1", "threshold"], ascending=[False, True]).iloc[0].threshold)\n', 'threshold_scores.to_csv(OUTPUT_ROOT / "roberta_validation_threshold_search.csv", index=False)\n', '\n', 'idx_cal, idx_tune = train_test_split(np.arange(len(val)), test_size=0.5, random_state=SEED, stratify=val.label)\n', 'def logit(p):\n', '    p = np.clip(np.asarray(p, float), 1e-6, 1-1e-6)\n', '    return np.log(p/(1-p)).reshape(-1,1)\n', 'platt = LogisticRegression(C=1e6, solver="lbfgs", random_state=SEED)\n', 'platt.fit(logit(val.p_text.iloc[idx_cal]), val.label.iloc[idx_cal])\n', 'p_tune = platt.predict_proba(logit(val.p_text.iloc[idx_tune]))[:,1]\n', 'platt_grid = pd.DataFrame({\n', '    "threshold": threshold_grid,\n', '    "tuning_half_macro_f1": [metrics(val.label.iloc[idx_tune], p_tune, t)["macro_f1"] for t in threshold_grid]\n', '})\n', 'platt_t = float(platt_grid.sort_values(["tuning_half_macro_f1", "threshold"], ascending=[False, True]).iloc[0].threshold)\n', 'platt_grid.to_csv(OUTPUT_ROOT / "roberta_platt_threshold_search.csv", index=False)\n', 'p_final_platt = platt.predict_proba(logit(final.probability_roberta))[:,1]\n', '\n', 'control_results = {\n', '    "roberta_default_0.5": metrics(final.label, final.probability_roberta, 0.5),\n', '    "roberta_validation_tuned_threshold": metrics(final.label, final.probability_roberta, best_t),\n', '    "roberta_platt_default_0.5": metrics(final.label, p_final_platt, 0.5),\n', '    "roberta_platt_tuned_threshold": metrics(final.label, p_final_platt, platt_t),\n', '    "locked_late_fusion": metrics(final.label, final.probability_fusion, 0.5),\n', '}\n', 'control_table = pd.DataFrame(control_results).T.reset_index(names="model")\n', 'control_table.to_csv(OUTPUT_ROOT / "fair_text_baseline_comparison.csv", index=False)\n', 'save_json("fair_text_baseline_comparison.json", {\n', '    "validation_selected_text_threshold": best_t,\n', '    "platt_calibration_fit_n": int(len(idx_cal)), "platt_threshold_tuning_n": int(len(idx_tune)),\n', '    "platt_selected_threshold": platt_t, "final_results": control_results\n', '})\n', 'display(control_table[["model","accuracy","macro_f1","roc_auc","pr_auc","brier","log_loss","threshold"]])']}, {'cell_type': 'markdown', 'id': '3ae0a2c3', 'metadata': {}, 'source': ['## 4. Source, domain, and time diagnostics\n', '\n', 'These are subgroup diagnostics, not a source-disjoint test: the trained models may have seen the same source categories during training. A source-only baseline is also fitted from original training labels. If it performs well, source identity alone carries target information and remains a plausible shortcut even though metadata was withheld from the neural networks.']}, {'cell_type': 'code', 'execution_count': None, 'id': '3d920cb2', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:58.611082Z', 'iopub.status.busy': '2026-09-09T12:46:58.611082Z', 'iopub.status.idle': '2026-09-09T12:47:00.701071Z', 'shell.execute_reply': '2026-09-09T12:47:00.701071Z'}}, 'outputs': [], 'source': ['test_meta = read_raw("test", ["id","subreddit","domain","created_utc","2_way_label"])\n', 'test_meta["id"] = test_meta["id"].astype(str); final["id"] = final["id"].astype(str)\n', 'enriched = final.merge(test_meta, on="id", how="left", validate="one_to_one")\n', 'enriched["year"] = pd.to_datetime(enriched.created_utc, unit="s", errors="coerce", utc=True).dt.year\n', '\n', 'def subgroup_table(group, min_n=30):\n', '    rows=[]\n', '    for key, g in enriched.groupby(group, dropna=False):\n', '        if len(g) < min_n or g.label.nunique() < 2: continue\n', '        tm=metrics(g.label, g.probability_roberta); fm=metrics(g.label, g.probability_fusion)\n', '        rows.append({group:key, "n":len(g), "class_1_rate":g.label.mean(),\n', '                     "roberta_macro_f1":tm["macro_f1"], "fusion_macro_f1":fm["macro_f1"],\n', '                     "fusion_delta_macro_f1":fm["macro_f1"]-tm["macro_f1"],\n', '                     "roberta_accuracy":tm["accuracy"], "fusion_accuracy":fm["accuracy"]})\n', '    columns=[group,"n","class_1_rate","roberta_macro_f1","fusion_macro_f1",\n', '             "fusion_delta_macro_f1","roberta_accuracy","fusion_accuracy"]\n', '    return pd.DataFrame(rows, columns=columns).sort_values("n", ascending=False)\n', '\n', 'for group in ["subreddit","domain","year"]:\n', '    table=subgroup_table(group)\n', '    table.to_csv(OUTPUT_ROOT / f"final_performance_by_{group}.csv", index=False)\n', '    display(table.head(15))\n', '\n', 'train_source = read_raw("train", ["subreddit","2_way_label"])\n', 'global_rate = float(train_source["2_way_label"].mean())\n', 'rates = train_source.groupby("subreddit")["2_way_label"].agg(["mean","size"])\n', 'smooth = (rates["mean"]*rates["size"] + global_rate*50)/(rates["size"]+50)\n', 'source_prob = enriched["subreddit"].map(smooth).fillna(global_rate).to_numpy()\n', 'source_only = metrics(enriched.label, source_prob, 0.5)\n', '\n', 'source_label_tab = pd.crosstab(train_source.subreddit, train_source["2_way_label"])\n', 'chi2, p, _, _ = chi2_contingency(source_label_tab)\n', 'v = math.sqrt(chi2/(source_label_tab.to_numpy().sum()*min(source_label_tab.shape[0]-1, source_label_tab.shape[1]-1)))\n', 'source_summary={"source_only_final_holdout":source_only,"training_source_label_cramers_v":float(v),"chi_square_p":float(p)}\n', 'save_json("source_shortcut_audit.json", source_summary)\n', 'print(source_summary)']}, {'cell_type': 'markdown', 'id': 'e1ded58e', 'metadata': {}, 'source': ['## 5. Perceptual duplicate screening\n', '\n', 'Exact hashes miss resized or recompressed copies. A 64-bit perceptual hash is computed for every usable development image and final image. A BK-tree searches for cross-set pairs within Hamming distance 6. These pairs are candidates for manual review; perceptual similarity alone is not proof of duplication.']}, {'cell_type': 'code', 'execution_count': None, 'id': '4ad4e1df', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:47:00.703077Z', 'iopub.status.busy': '2026-09-09T12:47:00.703077Z', 'iopub.status.idle': '2026-09-09T12:47:20.723448Z', 'shell.execute_reply': '2026-09-09T12:47:20.722944Z'}}, 'outputs': [], 'source': ['def resolve_original(path_value):\n', '    p=Path(str(path_value)); return p if p.is_absolute() else ORIGINAL_ROOT/p\n', '\n', 'def phash64(path):\n', '    with Image.open(path) as im:\n', '        a=np.asarray(im.convert("L").resize((32,32), Image.Resampling.LANCZOS), dtype=float)\n', '    low=dctn(a, type=2, norm="ortho")[:8,:8]\n', '    med=np.median(low.ravel()[1:])\n', '    bits=(low>med).ravel()\n', '    value=0\n', '    for bit in bits: value=(value<<1)|int(bit)\n', '    return value\n', '\n', 'cache_path=OUTPUT_ROOT/"perceptual_hashes.csv"\n', 'if cache_path.exists():\n', '    hashes=pd.read_csv(cache_path, dtype={"id":str,"phash_hex":str})\n', 'else:\n', '    image_rows=[]\n', '    for split in ["train","validation","test"]:\n', '        d=pd.read_parquet(PROCESSED_ROOT/"development_clean"/f"{split}.parquet")\n', '        image_rows.extend(("development",str(r.id),resolve_original(r.image_path)) for r in d.itertuples())\n', '    hold=pd.read_parquet(PROCESSED_ROOT/"final_holdout"/"final_5000.parquet")\n', '    image_rows.extend(("final",str(r.id),resolve_original(r.image_path)) for r in hold.itertuples())\n', '    out=[]\n', '    for i,(partition,sid,path) in enumerate(image_rows,1):\n', '        try: out.append({"partition":partition,"id":sid,"path":str(path),"phash_hex":f"{phash64(path):016x}","error":""})\n', '        except Exception as e: out.append({"partition":partition,"id":sid,"path":str(path),"phash_hex":"","error":type(e).__name__})\n', '        if i%2500==0: print(f"Hashed {i:,}/{len(image_rows):,}")\n', '    hashes=pd.DataFrame(out); hashes.to_csv(cache_path,index=False)\n', '\n', 'class BKNode:\n', '    def __init__(self,key,payload): self.key,self.payload,self.children=key,[payload],{}\n', '    def add(self,key,payload):\n', '        node=self\n', '        while True:\n', '            dist=(node.key^key).bit_count()\n', '            if dist==0: node.payload.append(payload); return\n', '            if dist not in node.children: node.children[dist]=BKNode(key,payload); return\n', '            node=node.children[dist]\n', '    def search(self,key,radius):\n', '        found=[]; stack=[self]\n', '        while stack:\n', '            node=stack.pop(); dist=(node.key^key).bit_count()\n', '            if dist<=radius: found.extend((p,dist) for p in node.payload)\n', '            stack.extend(child for edge,child in node.children.items() if dist-radius<=edge<=dist+radius)\n', '        return found\n', '\n', 'dev=hashes[(hashes.partition=="development") & hashes.phash_hex.ne("")]\n', 'fin=hashes[(hashes.partition=="final") & hashes.phash_hex.ne("")]\n', 'tree=None\n', 'for r in dev.itertuples():\n', '    key=int(r.phash_hex,16)\n', '    if tree is None: tree=BKNode(key,(r.id,r.path,r.phash_hex))\n', '    else: tree.add(key,(r.id,r.path,r.phash_hex))\n', 'pairs=[]\n', 'for r in fin.itertuples():\n', '    for (dev_id,dev_path,dev_hash),distance in tree.search(int(r.phash_hex,16),6):\n', '        pairs.append({"final_id":r.id,"development_id":dev_id,"hamming_distance":distance,\n', '                      "final_path":r.path,"development_path":dev_path,"final_phash":r.phash_hex,"development_phash":dev_hash})\n', 'near=pd.DataFrame(pairs).sort_values(["hamming_distance","final_id"]) if pairs else pd.DataFrame(columns=["final_id","development_id","hamming_distance"])\n', 'near.to_csv(OUTPUT_ROOT/"perceptual_near_duplicate_candidates.csv",index=False)\n', 'print(f"Usable hashes: development={len(dev):,}; final={len(fin):,}")\n', 'print(f"Cross-set candidate pairs at Hamming distance <=6: {len(near):,}")\n', 'display(near.head(20))']}, {'cell_type': 'markdown', 'id': 'ec90d45b', 'metadata': {}, 'source': ['## 6. Stronger split manifests for future retraining\n', '\n', 'The current checkpoints cannot be converted into source-disjoint or chronological experiments after training. This section creates reproducible manifests for those experiments without running expensive model training. Each manifest uses only the existing cleaned multimodal development examples.']}, {'cell_type': 'code', 'execution_count': None, 'id': '5a6267a2', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:47:20.726453Z', 'iopub.status.busy': '2026-09-09T12:47:20.725454Z', 'iopub.status.idle': '2026-09-09T12:47:24.549646Z', 'shell.execute_reply': '2026-09-09T12:47:24.549646Z'}}, 'outputs': [], 'source': ['clean_parts=[]\n', 'for split in ["train","validation","test"]:\n', '    d=pd.read_parquet(PROCESSED_ROOT/"development_clean"/f"{split}.parquet")\n', '    meta=read_raw(split,["id","subreddit","domain","created_utc","2_way_label"])\n', '    d["id"]=d.id.astype(str); meta["id"]=meta.id.astype(str)\n', '    clean_parts.append(d.merge(meta,on="id",how="left",validate="one_to_one"))\n', 'clean=pd.concat(clean_parts,ignore_index=True).drop_duplicates("id")\n', 'clean["created_datetime"]=pd.to_datetime(clean.created_utc,unit="s",errors="coerce",utc=True)\n', '\n', '# Source-disjoint: Fakeddit subreddits are label-pure. Allocate whole subreddits\n', '# separately inside each label so every split contains both classes.\n', 'purity=clean.groupby("subreddit")["label"].nunique()\n', 'assert purity.max()==1, "Expected subreddit-level distant-supervision labels."\n', 'source_labels=clean.groupby("subreddit")["label"].first()\n', 'counts=clean.groupby("subreddit").size()\n', 'assignment={}\n', 'for label in sorted(clean.label.unique()):\n', '    label_counts=counts[source_labels==label].sort_values(ascending=False)\n', '    label_total=int(label_counts.sum())\n', '    targets={"train":.70*label_total,"validation":.15*label_total,"test":.15*label_total}\n', '    totals={k:0 for k in targets}\n', '    for source,count in label_counts.items():\n', '        split=min(targets,key=lambda k: totals[k]/targets[k])\n', '        assignment[source]=split; totals[split]+=int(count)\n', 'source_manifest=clean[["id","label","text","image_path","subreddit","domain","created_utc"]].copy()\n', 'source_manifest["v2_split"]=source_manifest.subreddit.map(assignment)\n', 'assert source_manifest.groupby("subreddit").v2_split.nunique().max()==1\n', 'assert source_manifest.groupby("v2_split").label.nunique().min()==2\n', 'source_manifest.to_parquet(MANIFEST_ROOT/"source_disjoint.parquet",index=False)\n', '\n', 'chronological=clean.sort_values(["created_datetime","id"]).copy()\n', 'chronological["v2_split"]="train"\n', 'chronological.iloc[int(.70*len(chronological)):int(.85*len(chronological)), chronological.columns.get_loc("v2_split")]="validation"\n', 'chronological.iloc[int(.85*len(chronological)):, chronological.columns.get_loc("v2_split")]="test"\n', 'chronological[["id","label","text","image_path","subreddit","domain","created_utc","v2_split"]].to_parquet(\n', '    MANIFEST_ROOT/"chronological.parquet",index=False)\n', '\n', 'split_summary=pd.concat([\n', '    source_manifest.groupby("v2_split").agg(n=("id","size"),class_1_rate=("label","mean")).assign(manifest="source_disjoint"),\n', '    chronological.groupby("v2_split").agg(n=("id","size"),class_1_rate=("label","mean")).assign(manifest="chronological")\n', ']).reset_index()\n', 'split_summary.to_csv(OUTPUT_ROOT/"v2_manifest_summary.csv",index=False)\n', 'display(split_summary)']}, {'cell_type': 'markdown', 'id': '8d09aa3c', 'metadata': {}, 'source': ['## 7. Explainability coverage and reporting checks\n', '\n', 'This verifies whether the stored artifacts match the method description and writes a machine-readable correction list for the dissertation draft.']}, {'cell_type': 'code', 'execution_count': None, 'id': '9e0e1064', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:47:24.552126Z', 'iopub.status.busy': '2026-09-09T12:47:24.552126Z', 'iopub.status.idle': '2026-09-09T12:47:24.732109Z', 'shell.execute_reply': '2026-09-09T12:47:24.732109Z'}}, 'outputs': [], 'source': ['cases32=pd.read_csv(RESULTS_ROOT/"case_studies"/"all_32_multimodal_cases.csv")\n', 'cases8=pd.read_csv(RESULTS_ROOT/"case_studies"/"selected_8_case_studies.csv")\n', 'shap_summary=pd.read_csv(RESULTS_ROOT/"shap"/"shap_case_summary.csv")\n', 'grad_summary=pd.read_csv(RESULTS_ROOT/"gradcam"/"gradcam_case_summary.csv")\n', 'coverage={\n', '    "all_multimodal_cases":int(len(cases32)), "selected_paired_cases":int(len(cases8)),\n', '    "shap_cases":int(len(shap_summary)), "gradcam_cases":int(len(grad_summary)),\n', '    "case_columns":list(cases32.columns),\n', '}\n', 'if "label" in cases32.columns: coverage["all_32_label_counts"]={str(k):int(v) for k,v in cases32.label.value_counts().items()}\n', 'save_json("explainability_coverage.json",coverage)\n', '\n', 'raw_test_n=len(read_raw("test",["id"]))\n', 'robustness=json.loads((RESULTS_ROOT/"metrics"/"missing_modality_robustness"/"results.json").read_text())\n', 'changes={r["scenario"]:r["macro_f1_change_vs_full"] for r in robustness["results"]}\n', 'checks=pd.DataFrame([\n', '    {"item":"public test size","observed":raw_test_n,"expected":59319,"status":"PASS" if raw_test_n==59319 else "FAIL","draft_action":"Use 59,319 consistently."},\n', '    {"item":"missing text change sign","observed":changes.get("missing_text_image_fallback"),"expected":"negative","status":"PASS" if changes.get("missing_text_image_fallback",1)<0 else "FAIL","draft_action":"Report -0.0906, not +0.0906."},\n', '    {"item":"32-case table exists","observed":len(cases32),"expected":32,"status":"PASS" if len(cases32)==32 else "FAIL","draft_action":"Describe the full 32-case analysis and distinguish it from the four illustrated cases."},\n', '    {"item":"paired SHAP and Grad-CAM coverage","observed":f"SHAP={len(shap_summary)}, Grad-CAM={len(grad_summary)}","expected":">=32 each","status":"PASS" if min(len(shap_summary),len(grad_summary))>=32 else "FAIL","draft_action":"Reconcile claimed and generated explanation counts."},\n', '])\n', 'checks.to_csv(OUTPUT_ROOT/"reporting_consistency_checks.csv",index=False)\n', 'display(checks)\n', 'print(coverage)']}, {'cell_type': 'markdown', 'id': '2dda591b', 'metadata': {}, 'source': ['## Interpretation boundaries\n', '\n', 'The strongest supported conclusion remains specific: on the selected cleaned Fakeddit sample and locked checkpoints, late probability fusion improves over the original RoBERTa decision rule. The added controls show whether that advantage remains after fair threshold tuning and how strongly source and selection effects constrain generalisation.\n', '\n', 'The source-disjoint and chronological manifests must be used to retrain all models from scratch before making claims about transfer to unseen sources or later periods. Full training-seed uncertainty likewise requires several independent end-to-end training runs; it cannot be recovered from one checkpoint. This notebook deliberately does not fabricate those results.']}], 'metadata': {'kernelspec': {'display_name': 'Python 3', 'language': 'python', 'name': 'python3'}, 'language_info': {'codemirror_mode': {'name': 'ipython', 'version': 3}, 'file_extension': '.py', 'mimetype': 'text/x-python', 'name': 'python', 'nbconvert_exporter': 'python', 'pygments_lexer': 'ipython3', 'version': '3.12.3'}}, 'nbformat': 4, 'nbformat_minor': 5}, 'historical/v2/methodology_gap_analysis_v2.ipynb': {'cells': [{'cell_type': 'markdown', 'id': '4e390fca', 'metadata': {}, 'source': ['# Fakeddit multimodal methodology audit — v2\n', '\n', 'This notebook adds the methodological checks that were missing from the original project while preserving the original code, data, checkpoints, and results. It reads from `F:\\data sci\\project\\multimodal-fake-news-detection` and writes only to this `v2` folder.\n', '\n', 'The notebook covers:\n', '\n', '1. binary-label semantics and internal consistency;\n', '2. class-dependent image-selection bias;\n', '3. a fairer validation-tuned and calibrated RoBERTa comparison;\n', '4. source, domain, and time subgroup performance plus a source-only shortcut baseline;\n', '5. perceptual-image duplicate screening;\n', '6. source-disjoint and chronological manifests for stronger future retraining;\n', '7. explainability coverage and reporting consistency checks.\n', '\n', 'The final holdout is used only for locked evaluation of predeclared controls. No original model or result is overwritten.']}, {'cell_type': 'code', 'execution_count': 1, 'id': '150aecf6', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:48.042916Z', 'iopub.status.busy': '2026-09-09T12:46:48.041916Z', 'iopub.status.idle': '2026-09-09T12:46:49.845246Z', 'shell.execute_reply': '2026-09-09T12:46:49.845246Z'}}, 'outputs': [{'name': 'stdout', 'output_type': 'stream', 'text': ['Original (read-only): F:\\data sci\\project\\multimodal-fake-news-detection\n', 'v2 outputs: F:\\data sci\\project\\v2\n']}], 'source': ['from pathlib import Path\n', 'import json, hashlib, math, warnings\n', 'import numpy as np\n', 'import pandas as pd\n', 'import matplotlib.pyplot as plt\n', 'from PIL import Image\n', 'from scipy.fft import dctn\n', 'from scipy.stats import chi2_contingency\n', 'from sklearn.calibration import calibration_curve\n', 'from sklearn.linear_model import LogisticRegression\n', 'from sklearn.metrics import (\n', '    accuracy_score, precision_score, recall_score, f1_score,\n', '    roc_auc_score, average_precision_score, brier_score_loss,\n', '    log_loss, confusion_matrix\n', ')\n', 'from sklearn.model_selection import train_test_split\n', '\n', 'ORIGINAL_ROOT = Path(r"F:\\data sci\\project\\multimodal-fake-news-detection").resolve()\n', 'V2_ROOT = Path(r"F:\\data sci\\project\\v2").resolve()\n', 'OUTPUT_ROOT = V2_ROOT / "outputs"\n', 'MANIFEST_ROOT = V2_ROOT / "manifests"\n', 'RAW_ROOT = ORIGINAL_ROOT / "data" / "raw" / "fakeddit"\n', 'PROCESSED_ROOT = ORIGINAL_ROOT / "data" / "processed" / "fakeddit"\n', 'RESULTS_ROOT = ORIGINAL_ROOT / "results"\n', 'SEED = 2026\n', '\n', 'assert ORIGINAL_ROOT.exists(), ORIGINAL_ROOT\n', 'assert V2_ROOT != ORIGINAL_ROOT and ORIGINAL_ROOT not in V2_ROOT.parents\n', 'OUTPUT_ROOT.mkdir(parents=True, exist_ok=True)\n', 'MANIFEST_ROOT.mkdir(parents=True, exist_ok=True)\n', '\n', 'def save_json(name, obj):\n', '    path = OUTPUT_ROOT / name\n', '    path.write_text(json.dumps(obj, indent=2, default=str), encoding="utf-8")\n', '    return path\n', '\n', 'def raw_path(split):\n', '    name = {"train":"multimodal_train.tsv", "validation":"multimodal_validate.tsv", "test":"multimodal_test_public.tsv"}[split]\n', '    return RAW_ROOT / "multimodal_only_samples" / name\n', '\n', 'def read_raw(split, columns=None):\n', '    return pd.read_csv(raw_path(split), sep="\\t", usecols=columns, low_memory=False)\n', '\n', 'def metrics(y, p, threshold=0.5):\n', '    y = np.asarray(y, dtype=int); p = np.clip(np.asarray(p, dtype=float), 1e-7, 1-1e-7)\n', '    pred = (p >= threshold).astype(int)\n', '    return {\n', '        "n": int(len(y)), "threshold": float(threshold),\n', '        "accuracy": float(accuracy_score(y, pred)),\n', '        "precision": float(precision_score(y, pred, zero_division=0)),\n', '        "recall": float(recall_score(y, pred, zero_division=0)),\n', '        "f1": float(f1_score(y, pred, zero_division=0)),\n', '        "macro_f1": float(f1_score(y, pred, average="macro", zero_division=0)),\n', '        "roc_auc": float(roc_auc_score(y, p)) if len(np.unique(y)) == 2 else np.nan,\n', '        "pr_auc": float(average_precision_score(y, p)) if len(np.unique(y)) == 2 else np.nan,\n', '        "brier": float(brier_score_loss(y, p)),\n', '        "log_loss": float(log_loss(y, p, labels=[0,1])),\n', '        "confusion_matrix": confusion_matrix(y, pred, labels=[0,1]).tolist(),\n', '    }\n', '\n', 'print("Original (read-only):", ORIGINAL_ROOT)\n', 'print("v2 outputs:", V2_ROOT)']}, {'cell_type': 'markdown', 'id': '4d875460', 'metadata': {}, 'source': ['## 1. Verify label semantics\n', '\n', "Fakeddit's six-way label `0` is the true-content category; the other five categories are forms of false or misleading content. The binary encoding is therefore checked programmatically: binary class `1` must correspond exactly to six-way class `0`, and binary class `0` to six-way classes `1–5`."]}, {'cell_type': 'code', 'execution_count': 2, 'id': 'cf69b2b5', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:49.847787Z', 'iopub.status.busy': '2026-09-09T12:46:49.846782Z', 'iopub.status.idle': '2026-09-09T12:46:51.906215Z', 'shell.execute_reply': '2026-09-09T12:46:51.906215Z'}}, 'outputs': [{'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th>6_way_label</th>\n', '      <th>0</th>\n', '      <th>1</th>\n', '      <th>2</th>\n', '      <th>3</th>\n', '      <th>4</th>\n', '      <th>5</th>\n', '    </tr>\n', '    <tr>\n', '      <th>2_way_label</th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>0</td>\n', '      <td>33481</td>\n', '      <td>107221</td>\n', '      <td>11784</td>\n', '      <td>167857</td>\n', '      <td>21576</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>222081</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['6_way_label       0      1       2      3       4      5\n', '2_way_label                                             \n', '0                 0  33481  107221  11784  167857  21576\n', '1            222081      0       0      0       0      0']}, 'metadata': {}, 'output_type': 'display_data'}, {'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th>6_way_label</th>\n', '      <th>0</th>\n', '      <th>1</th>\n', '      <th>2</th>\n', '      <th>3</th>\n', '      <th>4</th>\n', '      <th>5</th>\n', '    </tr>\n', '    <tr>\n', '      <th>2_way_label</th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>0</td>\n', '      <td>3521</td>\n', '      <td>11277</td>\n', '      <td>1238</td>\n', '      <td>17810</td>\n', '      <td>2176</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>23320</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['6_way_label      0     1      2     3      4     5\n', '2_way_label                                       \n', '0                0  3521  11277  1238  17810  2176\n', '1            23320     0      0     0      0     0']}, 'metadata': {}, 'output_type': 'display_data'}, {'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th>6_way_label</th>\n', '      <th>0</th>\n', '      <th>1</th>\n', '      <th>2</th>\n', '      <th>3</th>\n', '      <th>4</th>\n', '      <th>5</th>\n', '    </tr>\n', '    <tr>\n', '      <th>2_way_label</th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '      <th></th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>0</td>\n', '      <td>3514</td>\n', '      <td>11297</td>\n', '      <td>1224</td>\n', '      <td>17472</td>\n', '      <td>2305</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>23507</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '      <td>0</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['6_way_label      0     1      2     3      4     5\n', '2_way_label                                       \n', '0                0  3514  11297  1224  17472  2305\n', '1            23507     0      0     0      0     0']}, 'metadata': {}, 'output_type': 'display_data'}, {'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>split</th>\n', '      <th>n</th>\n', '      <th>consistent_n</th>\n', '      <th>inconsistent_n</th>\n', '      <th>consistent_pct</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>train</td>\n', '      <td>564000</td>\n', '      <td>564000</td>\n', '      <td>0</td>\n', '      <td>100.0</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>validation</td>\n', '      <td>59342</td>\n', '      <td>59342</td>\n', '      <td>0</td>\n', '      <td>100.0</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>test</td>\n', '      <td>59319</td>\n', '      <td>59319</td>\n', '      <td>0</td>\n', '      <td>100.0</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['        split       n  consistent_n  inconsistent_n  consistent_pct\n', '0       train  564000        564000               0           100.0\n', '1  validation   59342         59342               0           100.0\n', '2        test   59319         59319               0           100.0']}, 'metadata': {}, 'output_type': 'display_data'}], 'source': ['label_rows = []\n', 'label_tables = {}\n', 'for split in ["train", "validation", "test"]:\n', '    d = read_raw(split, ["id", "2_way_label", "3_way_label", "6_way_label"])\n', '    tab = pd.crosstab(d["2_way_label"], d["6_way_label"])\n', '    label_tables[split] = tab\n', '    consistent = ((d["2_way_label"] == 1) == (d["6_way_label"] == 0))\n', '    label_rows.append({\n', '        "split": split, "n": len(d), "consistent_n": int(consistent.sum()),\n', '        "inconsistent_n": int((~consistent).sum()), "consistent_pct": float(100*consistent.mean())\n', '    })\n', '    display(tab)\n', '\n', 'label_audit = pd.DataFrame(label_rows)\n', 'label_audit.to_csv(OUTPUT_ROOT / "label_semantics_audit.csv", index=False)\n', 'assert label_audit["inconsistent_n"].sum() == 0\n', 'semantics = {\n', '    "binary_class_1": "true/real content",\n', '    "binary_class_0": "fake or misleading content (six-way classes 1-5)",\n', '    "verification": label_rows,\n', '    "limitation": "This verifies dataset encoding, not the factual correctness of every distant-supervision label."\n', '}\n', 'save_json("label_semantics.json", semantics)\n', 'display(label_audit)']}, {'cell_type': 'markdown', 'id': '3a8ba1ee', 'metadata': {}, 'source': ['## 2. Quantify selection bias caused by image availability\n', '\n', 'Equal sample IDs make comparisons between modalities fair within the retained subset. They do not make that subset representative. This section measures retention by label, year, domain, and subreddit and tests whether retention is independent of the binary label.']}, {'cell_type': 'code', 'execution_count': 3, 'id': 'de8fac17', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:51.908257Z', 'iopub.status.busy': '2026-09-09T12:46:51.908257Z', 'iopub.status.idle': '2026-09-09T12:46:55.460716Z', 'shell.execute_reply': '2026-09-09T12:46:55.460716Z'}}, 'outputs': [{'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>split</th>\n', '      <th>label</th>\n', '      <th>total</th>\n', '      <th>retained</th>\n', '      <th>retention_rate</th>\n', '      <th>removed</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>test</td>\n', '      <td>0</td>\n', '      <td>1811</td>\n', '      <td>861</td>\n', '      <td>0.475428</td>\n', '      <td>950</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>test</td>\n', '      <td>1</td>\n', '      <td>1189</td>\n', '      <td>1104</td>\n', '      <td>0.928511</td>\n', '      <td>85</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>train</td>\n', '      <td>0</td>\n', '      <td>12125</td>\n', '      <td>5854</td>\n', '      <td>0.482804</td>\n', '      <td>6271</td>\n', '    </tr>\n', '    <tr>\n', '      <th>3</th>\n', '      <td>train</td>\n', '      <td>1</td>\n', '      <td>7875</td>\n', '      <td>7275</td>\n', '      <td>0.923810</td>\n', '      <td>600</td>\n', '    </tr>\n', '    <tr>\n', '      <th>4</th>\n', '      <td>validation</td>\n', '      <td>0</td>\n', '      <td>1821</td>\n', '      <td>860</td>\n', '      <td>0.472268</td>\n', '      <td>961</td>\n', '    </tr>\n', '    <tr>\n', '      <th>5</th>\n', '      <td>validation</td>\n', '      <td>1</td>\n', '      <td>1179</td>\n', '      <td>1102</td>\n', '      <td>0.934690</td>\n', '      <td>77</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['        split  label  total  retained  retention_rate  removed\n', '0        test      0   1811       861        0.475428      950\n', '1        test      1   1189      1104        0.928511       85\n', '2       train      0  12125      5854        0.482804     6271\n', '3       train      1   7875      7275        0.923810      600\n', '4  validation      0   1821       860        0.472268      961\n', '5  validation      1   1179      1102        0.934690       77']}, 'metadata': {}, 'output_type': 'display_data'}, {'name': 'stdout', 'output_type': 'stream', 'text': ["{'n': 26000, 'chi_square': 5442.170120555753, 'p_value': 0.0, 'cramers_v': 0.4575087271364236, 'interpretation': 'Large dependence means complete-case filtering changes the target population. Macro-F1 does not remove this selection bias.'}\n"]}, {'data': {'image/png': '...', 'text/plain': ['<Figure size 700x400 with 1 Axes>']}, 'metadata': {}, 'output_type': 'display_data'}], 'source': ['status_parts = []\n', 'for split in ["train", "validation", "test"]:\n', '    p = PROCESSED_ROOT / "development_clean" / f"{split}_with_image_status.parquet"\n', '    s = pd.read_parquet(p)\n', '    meta = read_raw(split, ["id", "subreddit", "domain", "created_utc", "2_way_label"])\n', '    s["id"] = s["id"].astype(str); meta["id"] = meta["id"].astype(str)\n', '    s = s.merge(meta, on="id", how="left", validate="one_to_one")\n', '    s["retained"] = s["image_usable"].fillna(False).astype(bool)\n', '    s["year"] = pd.to_datetime(s["created_utc"], unit="s", errors="coerce", utc=True).dt.year\n', '    status_parts.append(s)\n', 'status = pd.concat(status_parts, ignore_index=True)\n', '\n', 'retention = (status.groupby(["split", "label"])["retained"]\n', '             .agg(total="size", retained="sum", retention_rate="mean").reset_index())\n', 'retention["removed"] = retention["total"] - retention["retained"]\n', 'retention.to_csv(OUTPUT_ROOT / "selection_retention_by_label.csv", index=False)\n', '\n', 'contingency = pd.crosstab(status["label"], status["retained"])\n', 'chi2, p_value, _, _ = chi2_contingency(contingency)\n', 'n = contingency.to_numpy().sum()\n', 'cramers_v = math.sqrt(chi2 / n)\n', 'bias_summary = {\n', '    "n": int(n), "chi_square": float(chi2), "p_value": float(p_value),\n', '    "cramers_v": float(cramers_v),\n', '    "interpretation": "Large dependence means complete-case filtering changes the target population. Macro-F1 does not remove this selection bias."\n', '}\n', 'save_json("selection_bias_summary.json", bias_summary)\n', '\n', 'for group in ["subreddit", "domain", "year"]:\n', '    g = (status.groupby(group, dropna=False)["retained"]\n', '         .agg(total="size", retained="sum", retention_rate="mean").reset_index())\n', '    g["removed"] = g["total"] - g["retained"]\n', '    g.sort_values(["total", "retention_rate"], ascending=[False, True]).to_csv(\n', '        OUTPUT_ROOT / f"selection_retention_by_{group}.csv", index=False)\n', '\n', 'display(retention)\n', 'print(bias_summary)\n', '\n', 'fig, ax = plt.subplots(figsize=(7,4))\n', 'for split, grp in retention.groupby("split"):\n', '    ax.plot(grp["label"].astype(str), grp["retention_rate"], marker="o", label=split)\n', 'ax.set(xlabel="Binary label (0=fake/misleading, 1=true)", ylabel="Image retention rate", ylim=(0,1),\n', '       title="Image filtering is strongly class-dependent")\n', 'ax.legend(); fig.tight_layout()\n', 'fig.savefig(OUTPUT_ROOT / "selection_retention_by_label.png", dpi=180)\n', 'plt.show()']}, {'cell_type': 'markdown', 'id': '0e54206c', 'metadata': {}, 'source': ['## 3. Fair text-only threshold and calibration controls\n', '\n', 'The original fusion weight was selected on validation macro-F1 while RoBERTa used the default 0.5 threshold. This section gives RoBERTa the same opportunity to tune its decision threshold. It also fits Platt calibration on one stratified half of validation and selects its threshold on the other half, then evaluates each predeclared variant once on the frozen holdout.']}, {'cell_type': 'code', 'execution_count': 4, 'id': '6fe2166a', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:55.462761Z', 'iopub.status.busy': '2026-09-09T12:46:55.462761Z', 'iopub.status.idle': '2026-09-09T12:46:58.608870Z', 'shell.execute_reply': '2026-09-09T12:46:58.608870Z'}}, 'outputs': [{'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>model</th>\n', '      <th>accuracy</th>\n', '      <th>macro_f1</th>\n', '      <th>roc_auc</th>\n', '      <th>pr_auc</th>\n', '      <th>brier</th>\n', '      <th>log_loss</th>\n', '      <th>threshold</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>roberta_default_0.5</td>\n', '      <td>0.8046</td>\n', '      <td>0.799966</td>\n', '      <td>0.884581</td>\n', '      <td>0.902735</td>\n', '      <td>0.151197</td>\n', '      <td>0.51234</td>\n', '      <td>0.5</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>roberta_validation_tuned_threshold</td>\n', '      <td>0.8038</td>\n', '      <td>0.800584</td>\n', '      <td>0.884581</td>\n', '      <td>0.902735</td>\n', '      <td>0.151197</td>\n', '      <td>0.51234</td>\n', '      <td>0.61</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>roberta_platt_default_0.5</td>\n', '      <td>0.805</td>\n', '      <td>0.800123</td>\n', '      <td>0.884581</td>\n', '      <td>0.902735</td>\n', '      <td>0.137634</td>\n', '      <td>0.430858</td>\n', '      <td>0.5</td>\n', '    </tr>\n', '    <tr>\n', '      <th>3</th>\n', '      <td>roberta_platt_tuned_threshold</td>\n', '      <td>0.8014</td>\n', '      <td>0.799667</td>\n', '      <td>0.884581</td>\n', '      <td>0.902735</td>\n', '      <td>0.137634</td>\n', '      <td>0.430858</td>\n', '      <td>0.64</td>\n', '    </tr>\n', '    <tr>\n', '      <th>4</th>\n', '      <td>locked_late_fusion</td>\n', '      <td>0.8242</td>\n', '      <td>0.818776</td>\n', '      <td>0.899306</td>\n', '      <td>0.909669</td>\n', '      <td>0.128115</td>\n', '      <td>0.404546</td>\n', '      <td>0.5</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['                                model accuracy  macro_f1   roc_auc    pr_auc  \\\n', '0                 roberta_default_0.5   0.8046  0.799966  0.884581  0.902735   \n', '1  roberta_validation_tuned_threshold   0.8038  0.800584  0.884581  0.902735   \n', '2           roberta_platt_default_0.5    0.805  0.800123  0.884581  0.902735   \n', '3       roberta_platt_tuned_threshold   0.8014  0.799667  0.884581  0.902735   \n', '4                  locked_late_fusion   0.8242  0.818776  0.899306  0.909669   \n', '\n', '      brier  log_loss threshold  \n', '0  0.151197   0.51234       0.5  \n', '1  0.151197   0.51234      0.61  \n', '2  0.137634  0.430858       0.5  \n', '3  0.137634  0.430858      0.64  \n', '4  0.128115  0.404546       0.5  ']}, 'metadata': {}, 'output_type': 'display_data'}], 'source': ['val = pd.read_csv(RESULTS_ROOT / "metrics" / "baseline_probabilities" / "roberta_validation.csv")\n', 'final = pd.read_csv(RESULTS_ROOT / "metrics" / "final_evaluation" / "final_predictions.csv")\n', 'val = val.rename(columns={"probability_class_1":"p_text"})\n', '\n', 'threshold_grid = np.linspace(0.05, 0.95, 181)\n', 'threshold_scores = pd.DataFrame({\n', '    "threshold": threshold_grid,\n', '    "validation_macro_f1": [metrics(val.label, val.p_text, t)["macro_f1"] for t in threshold_grid]\n', '})\n', 'best_t = float(threshold_scores.sort_values(["validation_macro_f1", "threshold"], ascending=[False, True]).iloc[0].threshold)\n', 'threshold_scores.to_csv(OUTPUT_ROOT / "roberta_validation_threshold_search.csv", index=False)\n', '\n', 'idx_cal, idx_tune = train_test_split(np.arange(len(val)), test_size=0.5, random_state=SEED, stratify=val.label)\n', 'def logit(p):\n', '    p = np.clip(np.asarray(p, float), 1e-6, 1-1e-6)\n', '    return np.log(p/(1-p)).reshape(-1,1)\n', 'platt = LogisticRegression(C=1e6, solver="lbfgs", random_state=SEED)\n', 'platt.fit(logit(val.p_text.iloc[idx_cal]), val.label.iloc[idx_cal])\n', 'p_tune = platt.predict_proba(logit(val.p_text.iloc[idx_tune]))[:,1]\n', 'platt_grid = pd.DataFrame({\n', '    "threshold": threshold_grid,\n', '    "tuning_half_macro_f1": [metrics(val.label.iloc[idx_tune], p_tune, t)["macro_f1"] for t in threshold_grid]\n', '})\n', 'platt_t = float(platt_grid.sort_values(["tuning_half_macro_f1", "threshold"], ascending=[False, True]).iloc[0].threshold)\n', 'platt_grid.to_csv(OUTPUT_ROOT / "roberta_platt_threshold_search.csv", index=False)\n', 'p_final_platt = platt.predict_proba(logit(final.probability_roberta))[:,1]\n', '\n', 'control_results = {\n', '    "roberta_default_0.5": metrics(final.label, final.probability_roberta, 0.5),\n', '    "roberta_validation_tuned_threshold": metrics(final.label, final.probability_roberta, best_t),\n', '    "roberta_platt_default_0.5": metrics(final.label, p_final_platt, 0.5),\n', '    "roberta_platt_tuned_threshold": metrics(final.label, p_final_platt, platt_t),\n', '    "locked_late_fusion": metrics(final.label, final.probability_fusion, 0.5),\n', '}\n', 'control_table = pd.DataFrame(control_results).T.reset_index(names="model")\n', 'control_table.to_csv(OUTPUT_ROOT / "fair_text_baseline_comparison.csv", index=False)\n', 'save_json("fair_text_baseline_comparison.json", {\n', '    "validation_selected_text_threshold": best_t,\n', '    "platt_calibration_fit_n": int(len(idx_cal)), "platt_threshold_tuning_n": int(len(idx_tune)),\n', '    "platt_selected_threshold": platt_t, "final_results": control_results\n', '})\n', 'display(control_table[["model","accuracy","macro_f1","roc_auc","pr_auc","brier","log_loss","threshold"]])']}, {'cell_type': 'markdown', 'id': '3ae0a2c3', 'metadata': {}, 'source': ['## 4. Source, domain, and time diagnostics\n', '\n', 'These are subgroup diagnostics, not a source-disjoint test: the trained models may have seen the same source categories during training. A source-only baseline is also fitted from original training labels. If it performs well, source identity alone carries target information and remains a plausible shortcut even though metadata was withheld from the neural networks.']}, {'cell_type': 'code', 'execution_count': 5, 'id': '3d920cb2', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:46:58.611082Z', 'iopub.status.busy': '2026-09-09T12:46:58.611082Z', 'iopub.status.idle': '2026-09-09T12:47:00.701071Z', 'shell.execute_reply': '2026-09-09T12:47:00.701071Z'}}, 'outputs': [{'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>subreddit</th>\n', '      <th>n</th>\n', '      <th>class_1_rate</th>\n', '      <th>roberta_macro_f1</th>\n', '      <th>fusion_macro_f1</th>\n', '      <th>fusion_delta_macro_f1</th>\n', '      <th>roberta_accuracy</th>\n', '      <th>fusion_accuracy</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['Empty DataFrame\n', 'Columns: [subreddit, n, class_1_rate, roberta_macro_f1, fusion_macro_f1, fusion_delta_macro_f1, roberta_accuracy, fusion_accuracy]\n', 'Index: []']}, 'metadata': {}, 'output_type': 'display_data'}, {'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>domain</th>\n', '      <th>n</th>\n', '      <th>class_1_rate</th>\n', '      <th>roberta_macro_f1</th>\n', '      <th>fusion_macro_f1</th>\n', '      <th>fusion_delta_macro_f1</th>\n', '      <th>roberta_accuracy</th>\n', '      <th>fusion_accuracy</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>i.redd.it</td>\n', '      <td>2094</td>\n', '      <td>0.521968</td>\n', '      <td>0.817583</td>\n', '      <td>0.840956</td>\n', '      <td>0.023373</td>\n', '      <td>0.819007</td>\n', '      <td>0.842407</td>\n', '    </tr>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>i.imgur.com</td>\n', '      <td>967</td>\n', '      <td>0.535677</td>\n', '      <td>0.769624</td>\n', '      <td>0.819925</td>\n', '      <td>0.050301</td>\n', '      <td>0.770424</td>\n', '      <td>0.821096</td>\n', '    </tr>\n', '    <tr>\n', '      <th>3</th>\n', '      <td>imgur.com</td>\n', '      <td>391</td>\n', '      <td>0.248082</td>\n', '      <td>0.746168</td>\n', '      <td>0.769084</td>\n', '      <td>0.022916</td>\n', '      <td>0.790281</td>\n', '      <td>0.803069</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>i.reddituploads.com</td>\n', '      <td>52</td>\n', '      <td>0.461538</td>\n', '      <td>0.787755</td>\n', '      <td>0.787755</td>\n', '      <td>0.000000</td>\n', '      <td>0.788462</td>\n', '      <td>0.788462</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['                domain     n  class_1_rate  roberta_macro_f1  fusion_macro_f1  \\\n', '1            i.redd.it  2094      0.521968          0.817583         0.840956   \n', '0          i.imgur.com   967      0.535677          0.769624         0.819925   \n', '3            imgur.com   391      0.248082          0.746168         0.769084   \n', '2  i.reddituploads.com    52      0.461538          0.787755         0.787755   \n', '\n', '   fusion_delta_macro_f1  roberta_accuracy  fusion_accuracy  \n', '1               0.023373          0.819007         0.842407  \n', '0               0.050301          0.770424         0.821096  \n', '3               0.022916          0.790281         0.803069  \n', '2               0.000000          0.788462         0.788462  ']}, 'metadata': {}, 'output_type': 'display_data'}, {'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>year</th>\n', '      <th>n</th>\n', '      <th>class_1_rate</th>\n', '      <th>roberta_macro_f1</th>\n', '      <th>fusion_macro_f1</th>\n', '      <th>fusion_delta_macro_f1</th>\n', '      <th>roberta_accuracy</th>\n', '      <th>fusion_accuracy</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>7</th>\n', '      <td>2019</td>\n', '      <td>1632</td>\n', '      <td>0.689338</td>\n', '      <td>0.788266</td>\n', '      <td>0.817526</td>\n', '      <td>0.029261</td>\n', '      <td>0.816789</td>\n', '      <td>0.845588</td>\n', '    </tr>\n', '    <tr>\n', '      <th>6</th>\n', '      <td>2018</td>\n', '      <td>894</td>\n', '      <td>0.346756</td>\n', '      <td>0.800649</td>\n', '      <td>0.801694</td>\n', '      <td>0.001045</td>\n', '      <td>0.806488</td>\n', '      <td>0.806488</td>\n', '    </tr>\n', '    <tr>\n', '      <th>5</th>\n', '      <td>2017</td>\n', '      <td>803</td>\n', '      <td>0.412204</td>\n', '      <td>0.781150</td>\n', '      <td>0.795535</td>\n', '      <td>0.014385</td>\n', '      <td>0.782067</td>\n', '      <td>0.795766</td>\n', '    </tr>\n', '    <tr>\n', '      <th>4</th>\n', '      <td>2016</td>\n', '      <td>516</td>\n', '      <td>0.548450</td>\n', '      <td>0.805636</td>\n', '      <td>0.814241</td>\n', '      <td>0.008605</td>\n', '      <td>0.810078</td>\n', '      <td>0.819767</td>\n', '    </tr>\n', '    <tr>\n', '      <th>3</th>\n', '      <td>2015</td>\n', '      <td>434</td>\n', '      <td>0.640553</td>\n', '      <td>0.821607</td>\n', '      <td>0.821714</td>\n', '      <td>0.000107</td>\n', '      <td>0.836406</td>\n', '      <td>0.838710</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>2014</td>\n', '      <td>341</td>\n', '      <td>0.700880</td>\n', '      <td>0.739542</td>\n', '      <td>0.795830</td>\n', '      <td>0.056289</td>\n', '      <td>0.771261</td>\n', '      <td>0.821114</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>2013</td>\n', '      <td>240</td>\n', '      <td>0.633333</td>\n', '      <td>0.793681</td>\n', '      <td>0.836160</td>\n', '      <td>0.042478</td>\n', '      <td>0.800000</td>\n', '      <td>0.841667</td>\n', '    </tr>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>2012</td>\n', '      <td>127</td>\n', '      <td>0.606299</td>\n', '      <td>0.762587</td>\n', '      <td>0.801376</td>\n', '      <td>0.038789</td>\n', '      <td>0.763780</td>\n', '      <td>0.803150</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['   year     n  class_1_rate  roberta_macro_f1  fusion_macro_f1  \\\n', '7  2019  1632      0.689338          0.788266         0.817526   \n', '6  2018   894      0.346756          0.800649         0.801694   \n', '5  2017   803      0.412204          0.781150         0.795535   \n', '4  2016   516      0.548450          0.805636         0.814241   \n', '3  2015   434      0.640553          0.821607         0.821714   \n', '2  2014   341      0.700880          0.739542         0.795830   \n', '1  2013   240      0.633333          0.793681         0.836160   \n', '0  2012   127      0.606299          0.762587         0.801376   \n', '\n', '   fusion_delta_macro_f1  roberta_accuracy  fusion_accuracy  \n', '7               0.029261          0.816789         0.845588  \n', '6               0.001045          0.806488         0.806488  \n', '5               0.014385          0.782067         0.795766  \n', '4               0.008605          0.810078         0.819767  \n', '3               0.000107          0.836406         0.838710  \n', '2               0.056289          0.771261         0.821114  \n', '1               0.042478          0.800000         0.841667  \n', '0               0.038789          0.763780         0.803150  ']}, 'metadata': {}, 'output_type': 'display_data'}, {'name': 'stdout', 'output_type': 'stream', 'text': ["{'source_only_final_holdout': {'n': 5000, 'threshold': 0.5, 'accuracy': 1.0, 'precision': 1.0, 'recall': 1.0, 'f1': 1.0, 'macro_f1': 1.0, 'roc_auc': 0.9999999999999999, 'pr_auc': 1.0, 'brier': 8.307496693354844e-06, 'log_loss': 0.0012454003788193238, 'confusion_matrix': [[2201, 0], [0, 2799]]}, 'training_source_label_cramers_v': 1.0, 'chi_square_p': 0.0}\n"]}], 'source': ['test_meta = read_raw("test", ["id","subreddit","domain","created_utc","2_way_label"])\n', 'test_meta["id"] = test_meta["id"].astype(str); final["id"] = final["id"].astype(str)\n', 'enriched = final.merge(test_meta, on="id", how="left", validate="one_to_one")\n', 'enriched["year"] = pd.to_datetime(enriched.created_utc, unit="s", errors="coerce", utc=True).dt.year\n', '\n', 'def subgroup_table(group, min_n=30):\n', '    rows=[]\n', '    for key, g in enriched.groupby(group, dropna=False):\n', '        if len(g) < min_n or g.label.nunique() < 2: continue\n', '        tm=metrics(g.label, g.probability_roberta); fm=metrics(g.label, g.probability_fusion)\n', '        rows.append({group:key, "n":len(g), "class_1_rate":g.label.mean(),\n', '                     "roberta_macro_f1":tm["macro_f1"], "fusion_macro_f1":fm["macro_f1"],\n', '                     "fusion_delta_macro_f1":fm["macro_f1"]-tm["macro_f1"],\n', '                     "roberta_accuracy":tm["accuracy"], "fusion_accuracy":fm["accuracy"]})\n', '    columns=[group,"n","class_1_rate","roberta_macro_f1","fusion_macro_f1",\n', '             "fusion_delta_macro_f1","roberta_accuracy","fusion_accuracy"]\n', '    return pd.DataFrame(rows, columns=columns).sort_values("n", ascending=False)\n', '\n', 'for group in ["subreddit","domain","year"]:\n', '    table=subgroup_table(group)\n', '    table.to_csv(OUTPUT_ROOT / f"final_performance_by_{group}.csv", index=False)\n', '    display(table.head(15))\n', '\n', 'train_source = read_raw("train", ["subreddit","2_way_label"])\n', 'global_rate = float(train_source["2_way_label"].mean())\n', 'rates = train_source.groupby("subreddit")["2_way_label"].agg(["mean","size"])\n', 'smooth = (rates["mean"]*rates["size"] + global_rate*50)/(rates["size"]+50)\n', 'source_prob = enriched["subreddit"].map(smooth).fillna(global_rate).to_numpy()\n', 'source_only = metrics(enriched.label, source_prob, 0.5)\n', '\n', 'source_label_tab = pd.crosstab(train_source.subreddit, train_source["2_way_label"])\n', 'chi2, p, _, _ = chi2_contingency(source_label_tab)\n', 'v = math.sqrt(chi2/(source_label_tab.to_numpy().sum()*min(source_label_tab.shape[0]-1, source_label_tab.shape[1]-1)))\n', 'source_summary={"source_only_final_holdout":source_only,"training_source_label_cramers_v":float(v),"chi_square_p":float(p)}\n', 'save_json("source_shortcut_audit.json", source_summary)\n', 'print(source_summary)']}, {'cell_type': 'markdown', 'id': 'e1ded58e', 'metadata': {}, 'source': ['## 5. Perceptual duplicate screening\n', '\n', 'Exact hashes miss resized or recompressed copies. A 64-bit perceptual hash is computed for every usable development image and final image. A BK-tree searches for cross-set pairs within Hamming distance 6. These pairs are candidates for manual review; perceptual similarity alone is not proof of duplication.']}, {'cell_type': 'code', 'execution_count': 6, 'id': '4ad4e1df', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:47:00.703077Z', 'iopub.status.busy': '2026-09-09T12:47:00.703077Z', 'iopub.status.idle': '2026-09-09T12:47:20.723448Z', 'shell.execute_reply': '2026-09-09T12:47:20.722944Z'}}, 'outputs': [{'name': 'stdout', 'output_type': 'stream', 'text': ['Usable hashes: development=17,056; final=5,000\n', 'Cross-set candidate pairs at Hamming distance <=6: 45\n']}, {'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>final_id</th>\n', '      <th>development_id</th>\n', '      <th>hamming_distance</th>\n', '      <th>final_path</th>\n', '      <th>development_path</th>\n', '      <th>final_phash</th>\n', '      <th>development_phash</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>36</th>\n', '      <td>1f7ss5</td>\n', '      <td>22gc0g</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>87c330e535da6b0d</td>\n', '      <td>87c330e535da6b0d</td>\n', '    </tr>\n', '    <tr>\n', '      <th>13</th>\n', '      <td>1nyf1b</td>\n', '      <td>1nv0il</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>ee4743131e3e36a1</td>\n', '      <td>ee4743131e3e36a1</td>\n', '    </tr>\n', '    <tr>\n', '      <th>10</th>\n', '      <td>1utjen</td>\n', '      <td>5q44vv</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>d2342fca70c3ce9c</td>\n', '      <td>d2342fca70c3ce9c</td>\n', '    </tr>\n', '    <tr>\n', '      <th>11</th>\n', '      <td>1utjen</td>\n', '      <td>5z7g98</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>d2342fca70c3ce9c</td>\n', '      <td>d2342fca70c3ce9c</td>\n', '    </tr>\n', '    <tr>\n', '      <th>12</th>\n', '      <td>1utjen</td>\n', '      <td>3gzmch</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>d2342fca70c3ce9c</td>\n', '      <td>d2342fca70c3ce9c</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>2mzoha</td>\n', '      <td>azf49b</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>efc5903ab2644d8d</td>\n', '      <td>efc5903ab2644d8d</td>\n', '    </tr>\n', '    <tr>\n', '      <th>32</th>\n', '      <td>3pi4te</td>\n', '      <td>5wpg4c</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>9209ab3e3cd86aa7</td>\n', '      <td>9209ab3e3cd86aa7</td>\n', '    </tr>\n', '    <tr>\n', '      <th>19</th>\n', '      <td>4naxwc</td>\n', '      <td>51qjm4</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>8000000000000000</td>\n', '      <td>8000000000000000</td>\n', '    </tr>\n', '    <tr>\n', '      <th>20</th>\n', '      <td>4naxwc</td>\n', '      <td>7uv14s</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>8000000000000000</td>\n', '      <td>8000000000000000</td>\n', '    </tr>\n', '    <tr>\n', '      <th>21</th>\n', '      <td>4naxwc</td>\n', '      <td>cw2u0g</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>8000000000000000</td>\n', '      <td>8000000000000000</td>\n', '    </tr>\n', '    <tr>\n', '      <th>22</th>\n', '      <td>4naxwc</td>\n', '      <td>chab3g</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>8000000000000000</td>\n', '      <td>8000000000000000</td>\n', '    </tr>\n', '    <tr>\n', '      <th>23</th>\n', '      <td>4naxwc</td>\n', '      <td>cyt4eo</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>8000000000000000</td>\n', '      <td>8000000000000000</td>\n', '    </tr>\n', '    <tr>\n', '      <th>24</th>\n', '      <td>4naxwc</td>\n', '      <td>8my9h0</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>8000000000000000</td>\n', '      <td>8000000000000000</td>\n', '    </tr>\n', '    <tr>\n', '      <th>14</th>\n', '      <td>4snxdo</td>\n', '      <td>25dl0y</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>b682f2309e26e71e</td>\n', '      <td>b682f2309e26e71e</td>\n', '    </tr>\n', '    <tr>\n', '      <th>42</th>\n', '      <td>4wwwx1</td>\n', '      <td>4icuhx</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>c0c0c060ecfeeef9</td>\n', '      <td>c0c0c060ecfeeef9</td>\n', '    </tr>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>50njnc</td>\n', '      <td>552nde</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>d03f2fd03b2fc0b0</td>\n', '      <td>d03f2fd03b2fc0b0</td>\n', '    </tr>\n', '    <tr>\n', '      <th>27</th>\n', '      <td>5htie8</td>\n', '      <td>75ccj4</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>f25a78b255f46289</td>\n', '      <td>f25a78b255f46289</td>\n', '    </tr>\n', '    <tr>\n', '      <th>44</th>\n', '      <td>6xep1b</td>\n', '      <td>9ewm59</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>d40f0fe7941f5813</td>\n', '      <td>d40f0fe7941f5813</td>\n', '    </tr>\n', '    <tr>\n', '      <th>26</th>\n', '      <td>7ce3a4</td>\n', '      <td>888xos</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>a06b5ada5a7c6616</td>\n', '      <td>a06b5ada5a7c6616</td>\n', '    </tr>\n', '    <tr>\n', '      <th>40</th>\n', '      <td>7frcnd</td>\n', '      <td>2zgjms</td>\n', '      <td>0</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>F:\\data sci\\project\\multimodal-fake-news-detec...</td>\n', '      <td>d44cec707237d613</td>\n', '      <td>d44cec707237d613</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['   final_id development_id  hamming_distance  \\\n', '36   1f7ss5         22gc0g                 0   \n', '13   1nyf1b         1nv0il                 0   \n', '10   1utjen         5q44vv                 0   \n', '11   1utjen         5z7g98                 0   \n', '12   1utjen         3gzmch                 0   \n', '1    2mzoha         azf49b                 0   \n', '32   3pi4te         5wpg4c                 0   \n', '19   4naxwc         51qjm4                 0   \n', '20   4naxwc         7uv14s                 0   \n', '21   4naxwc         cw2u0g                 0   \n', '22   4naxwc         chab3g                 0   \n', '23   4naxwc         cyt4eo                 0   \n', '24   4naxwc         8my9h0                 0   \n', '14   4snxdo         25dl0y                 0   \n', '42   4wwwx1         4icuhx                 0   \n', '0    50njnc         552nde                 0   \n', '27   5htie8         75ccj4                 0   \n', '44   6xep1b         9ewm59                 0   \n', '26   7ce3a4         888xos                 0   \n', '40   7frcnd         2zgjms                 0   \n', '\n', '                                           final_path  \\\n', '36  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '13  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '10  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '11  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '12  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '1   F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '32  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '19  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '20  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '21  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '22  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '23  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '24  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '14  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '42  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '0   F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '27  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '44  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '26  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '40  F:\\data sci\\project\\multimodal-fake-news-detec...   \n', '\n', '                                     development_path       final_phash  \\\n', '36  F:\\data sci\\project\\multimodal-fake-news-detec...  87c330e535da6b0d   \n', '13  F:\\data sci\\project\\multimodal-fake-news-detec...  ee4743131e3e36a1   \n', '10  F:\\data sci\\project\\multimodal-fake-news-detec...  d2342fca70c3ce9c   \n', '11  F:\\data sci\\project\\multimodal-fake-news-detec...  d2342fca70c3ce9c   \n', '12  F:\\data sci\\project\\multimodal-fake-news-detec...  d2342fca70c3ce9c   \n', '1   F:\\data sci\\project\\multimodal-fake-news-detec...  efc5903ab2644d8d   \n', '32  F:\\data sci\\project\\multimodal-fake-news-detec...  9209ab3e3cd86aa7   \n', '19  F:\\data sci\\project\\multimodal-fake-news-detec...  8000000000000000   \n', '20  F:\\data sci\\project\\multimodal-fake-news-detec...  8000000000000000   \n', '21  F:\\data sci\\project\\multimodal-fake-news-detec...  8000000000000000   \n', '22  F:\\data sci\\project\\multimodal-fake-news-detec...  8000000000000000   \n', '23  F:\\data sci\\project\\multimodal-fake-news-detec...  8000000000000000   \n', '24  F:\\data sci\\project\\multimodal-fake-news-detec...  8000000000000000   \n', '14  F:\\data sci\\project\\multimodal-fake-news-detec...  b682f2309e26e71e   \n', '42  F:\\data sci\\project\\multimodal-fake-news-detec...  c0c0c060ecfeeef9   \n', '0   F:\\data sci\\project\\multimodal-fake-news-detec...  d03f2fd03b2fc0b0   \n', '27  F:\\data sci\\project\\multimodal-fake-news-detec...  f25a78b255f46289   \n', '44  F:\\data sci\\project\\multimodal-fake-news-detec...  d40f0fe7941f5813   \n', '26  F:\\data sci\\project\\multimodal-fake-news-detec...  a06b5ada5a7c6616   \n', '40  F:\\data sci\\project\\multimodal-fake-news-detec...  d44cec707237d613   \n', '\n', '   development_phash  \n', '36  87c330e535da6b0d  \n', '13  ee4743131e3e36a1  \n', '10  d2342fca70c3ce9c  \n', '11  d2342fca70c3ce9c  \n', '12  d2342fca70c3ce9c  \n', '1   efc5903ab2644d8d  \n', '32  9209ab3e3cd86aa7  \n', '19  8000000000000000  \n', '20  8000000000000000  \n', '21  8000000000000000  \n', '22  8000000000000000  \n', '23  8000000000000000  \n', '24  8000000000000000  \n', '14  b682f2309e26e71e  \n', '42  c0c0c060ecfeeef9  \n', '0   d03f2fd03b2fc0b0  \n', '27  f25a78b255f46289  \n', '44  d40f0fe7941f5813  \n', '26  a06b5ada5a7c6616  \n', '40  d44cec707237d613  ']}, 'metadata': {}, 'output_type': 'display_data'}], 'source': ['def resolve_original(path_value):\n', '    p=Path(str(path_value)); return p if p.is_absolute() else ORIGINAL_ROOT/p\n', '\n', 'def phash64(path):\n', '    with Image.open(path) as im:\n', '        a=np.asarray(im.convert("L").resize((32,32), Image.Resampling.LANCZOS), dtype=float)\n', '    low=dctn(a, type=2, norm="ortho")[:8,:8]\n', '    med=np.median(low.ravel()[1:])\n', '    bits=(low>med).ravel()\n', '    value=0\n', '    for bit in bits: value=(value<<1)|int(bit)\n', '    return value\n', '\n', 'cache_path=OUTPUT_ROOT/"perceptual_hashes.csv"\n', 'if cache_path.exists():\n', '    hashes=pd.read_csv(cache_path, dtype={"id":str,"phash_hex":str})\n', 'else:\n', '    image_rows=[]\n', '    for split in ["train","validation","test"]:\n', '        d=pd.read_parquet(PROCESSED_ROOT/"development_clean"/f"{split}.parquet")\n', '        image_rows.extend(("development",str(r.id),resolve_original(r.image_path)) for r in d.itertuples())\n', '    hold=pd.read_parquet(PROCESSED_ROOT/"final_holdout"/"final_5000.parquet")\n', '    image_rows.extend(("final",str(r.id),resolve_original(r.image_path)) for r in hold.itertuples())\n', '    out=[]\n', '    for i,(partition,sid,path) in enumerate(image_rows,1):\n', '        try: out.append({"partition":partition,"id":sid,"path":str(path),"phash_hex":f"{phash64(path):016x}","error":""})\n', '        except Exception as e: out.append({"partition":partition,"id":sid,"path":str(path),"phash_hex":"","error":type(e).__name__})\n', '        if i%2500==0: print(f"Hashed {i:,}/{len(image_rows):,}")\n', '    hashes=pd.DataFrame(out); hashes.to_csv(cache_path,index=False)\n', '\n', 'class BKNode:\n', '    def __init__(self,key,payload): self.key,self.payload,self.children=key,[payload],{}\n', '    def add(self,key,payload):\n', '        node=self\n', '        while True:\n', '            dist=(node.key^key).bit_count()\n', '            if dist==0: node.payload.append(payload); return\n', '            if dist not in node.children: node.children[dist]=BKNode(key,payload); return\n', '            node=node.children[dist]\n', '    def search(self,key,radius):\n', '        found=[]; stack=[self]\n', '        while stack:\n', '            node=stack.pop(); dist=(node.key^key).bit_count()\n', '            if dist<=radius: found.extend((p,dist) for p in node.payload)\n', '            stack.extend(child for edge,child in node.children.items() if dist-radius<=edge<=dist+radius)\n', '        return found\n', '\n', 'dev=hashes[(hashes.partition=="development") & hashes.phash_hex.ne("")]\n', 'fin=hashes[(hashes.partition=="final") & hashes.phash_hex.ne("")]\n', 'tree=None\n', 'for r in dev.itertuples():\n', '    key=int(r.phash_hex,16)\n', '    if tree is None: tree=BKNode(key,(r.id,r.path,r.phash_hex))\n', '    else: tree.add(key,(r.id,r.path,r.phash_hex))\n', 'pairs=[]\n', 'for r in fin.itertuples():\n', '    for (dev_id,dev_path,dev_hash),distance in tree.search(int(r.phash_hex,16),6):\n', '        pairs.append({"final_id":r.id,"development_id":dev_id,"hamming_distance":distance,\n', '                      "final_path":r.path,"development_path":dev_path,"final_phash":r.phash_hex,"development_phash":dev_hash})\n', 'near=pd.DataFrame(pairs).sort_values(["hamming_distance","final_id"]) if pairs else pd.DataFrame(columns=["final_id","development_id","hamming_distance"])\n', 'near.to_csv(OUTPUT_ROOT/"perceptual_near_duplicate_candidates.csv",index=False)\n', 'print(f"Usable hashes: development={len(dev):,}; final={len(fin):,}")\n', 'print(f"Cross-set candidate pairs at Hamming distance <=6: {len(near):,}")\n', 'display(near.head(20))']}, {'cell_type': 'markdown', 'id': 'ec90d45b', 'metadata': {}, 'source': ['## 6. Stronger split manifests for future retraining\n', '\n', 'The current checkpoints cannot be converted into source-disjoint or chronological experiments after training. This section creates reproducible manifests for those experiments without running expensive model training. Each manifest uses only the existing cleaned multimodal development examples.']}, {'cell_type': 'code', 'execution_count': 7, 'id': '5a6267a2', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:47:20.726453Z', 'iopub.status.busy': '2026-09-09T12:47:20.725454Z', 'iopub.status.idle': '2026-09-09T12:47:24.549646Z', 'shell.execute_reply': '2026-09-09T12:47:24.549646Z'}}, 'outputs': [{'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>v2_split</th>\n', '      <th>n</th>\n', '      <th>class_1_rate</th>\n', '      <th>manifest</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>test</td>\n', '      <td>2739</td>\n', '      <td>0.546915</td>\n', '      <td>source_disjoint</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>train</td>\n', '      <td>10524</td>\n', '      <td>0.529171</td>\n', '      <td>source_disjoint</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>validation</td>\n', '      <td>3793</td>\n', '      <td>0.636436</td>\n', '      <td>source_disjoint</td>\n', '    </tr>\n', '    <tr>\n', '      <th>3</th>\n', '      <td>test</td>\n', '      <td>2559</td>\n', '      <td>0.711606</td>\n', '      <td>chronological</td>\n', '    </tr>\n', '    <tr>\n', '      <th>4</th>\n', '      <td>train</td>\n', '      <td>11939</td>\n', '      <td>0.500377</td>\n', '      <td>chronological</td>\n', '    </tr>\n', '    <tr>\n', '      <th>5</th>\n', '      <td>validation</td>\n', '      <td>2558</td>\n', '      <td>0.659109</td>\n', '      <td>chronological</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['     v2_split      n  class_1_rate         manifest\n', '0        test   2739      0.546915  source_disjoint\n', '1       train  10524      0.529171  source_disjoint\n', '2  validation   3793      0.636436  source_disjoint\n', '3        test   2559      0.711606    chronological\n', '4       train  11939      0.500377    chronological\n', '5  validation   2558      0.659109    chronological']}, 'metadata': {}, 'output_type': 'display_data'}], 'source': ['clean_parts=[]\n', 'for split in ["train","validation","test"]:\n', '    d=pd.read_parquet(PROCESSED_ROOT/"development_clean"/f"{split}.parquet")\n', '    meta=read_raw(split,["id","subreddit","domain","created_utc","2_way_label"])\n', '    d["id"]=d.id.astype(str); meta["id"]=meta.id.astype(str)\n', '    clean_parts.append(d.merge(meta,on="id",how="left",validate="one_to_one"))\n', 'clean=pd.concat(clean_parts,ignore_index=True).drop_duplicates("id")\n', 'clean["created_datetime"]=pd.to_datetime(clean.created_utc,unit="s",errors="coerce",utc=True)\n', '\n', '# Source-disjoint: Fakeddit subreddits are label-pure. Allocate whole subreddits\n', '# separately inside each label so every split contains both classes.\n', 'purity=clean.groupby("subreddit")["label"].nunique()\n', 'assert purity.max()==1, "Expected subreddit-level distant-supervision labels."\n', 'source_labels=clean.groupby("subreddit")["label"].first()\n', 'counts=clean.groupby("subreddit").size()\n', 'assignment={}\n', 'for label in sorted(clean.label.unique()):\n', '    label_counts=counts[source_labels==label].sort_values(ascending=False)\n', '    label_total=int(label_counts.sum())\n', '    targets={"train":.70*label_total,"validation":.15*label_total,"test":.15*label_total}\n', '    totals={k:0 for k in targets}\n', '    for source,count in label_counts.items():\n', '        split=min(targets,key=lambda k: totals[k]/targets[k])\n', '        assignment[source]=split; totals[split]+=int(count)\n', 'source_manifest=clean[["id","label","text","image_path","subreddit","domain","created_utc"]].copy()\n', 'source_manifest["v2_split"]=source_manifest.subreddit.map(assignment)\n', 'assert source_manifest.groupby("subreddit").v2_split.nunique().max()==1\n', 'assert source_manifest.groupby("v2_split").label.nunique().min()==2\n', 'source_manifest.to_parquet(MANIFEST_ROOT/"source_disjoint.parquet",index=False)\n', '\n', 'chronological=clean.sort_values(["created_datetime","id"]).copy()\n', 'chronological["v2_split"]="train"\n', 'chronological.iloc[int(.70*len(chronological)):int(.85*len(chronological)), chronological.columns.get_loc("v2_split")]="validation"\n', 'chronological.iloc[int(.85*len(chronological)):, chronological.columns.get_loc("v2_split")]="test"\n', 'chronological[["id","label","text","image_path","subreddit","domain","created_utc","v2_split"]].to_parquet(\n', '    MANIFEST_ROOT/"chronological.parquet",index=False)\n', '\n', 'split_summary=pd.concat([\n', '    source_manifest.groupby("v2_split").agg(n=("id","size"),class_1_rate=("label","mean")).assign(manifest="source_disjoint"),\n', '    chronological.groupby("v2_split").agg(n=("id","size"),class_1_rate=("label","mean")).assign(manifest="chronological")\n', ']).reset_index()\n', 'split_summary.to_csv(OUTPUT_ROOT/"v2_manifest_summary.csv",index=False)\n', 'display(split_summary)']}, {'cell_type': 'markdown', 'id': '8d09aa3c', 'metadata': {}, 'source': ['## 7. Explainability coverage and reporting checks\n', '\n', 'This verifies whether the stored artifacts match the method description and writes a machine-readable correction list for the dissertation draft.']}, {'cell_type': 'code', 'execution_count': 8, 'id': '9e0e1064', 'metadata': {'execution': {'iopub.execute_input': '2026-09-09T12:47:24.552126Z', 'iopub.status.busy': '2026-09-09T12:47:24.552126Z', 'iopub.status.idle': '2026-09-09T12:47:24.732109Z', 'shell.execute_reply': '2026-09-09T12:47:24.732109Z'}}, 'outputs': [{'data': {'text/html': ['<div>\n', '<style scoped>\n', '    .dataframe tbody tr th:only-of-type {\n', '        vertical-align: middle;\n', '    }\n', '\n', '    .dataframe tbody tr th {\n', '        vertical-align: top;\n', '    }\n', '\n', '    .dataframe thead th {\n', '        text-align: right;\n', '    }\n', '</style>\n', '<table border="1" class="dataframe">\n', '  <thead>\n', '    <tr style="text-align: right;">\n', '      <th></th>\n', '      <th>item</th>\n', '      <th>observed</th>\n', '      <th>expected</th>\n', '      <th>status</th>\n', '      <th>draft_action</th>\n', '    </tr>\n', '  </thead>\n', '  <tbody>\n', '    <tr>\n', '      <th>0</th>\n', '      <td>public test size</td>\n', '      <td>59319</td>\n', '      <td>59319</td>\n', '      <td>PASS</td>\n', '      <td>Use 59,319 consistently.</td>\n', '    </tr>\n', '    <tr>\n', '      <th>1</th>\n', '      <td>missing text change sign</td>\n', '      <td>-0.090556</td>\n', '      <td>negative</td>\n', '      <td>PASS</td>\n', '      <td>Report -0.0906, not +0.0906.</td>\n', '    </tr>\n', '    <tr>\n', '      <th>2</th>\n', '      <td>32-case table exists</td>\n', '      <td>32</td>\n', '      <td>32</td>\n', '      <td>PASS</td>\n', '      <td>Describe the full 32-case analysis and disting...</td>\n', '    </tr>\n', '    <tr>\n', '      <th>3</th>\n', '      <td>paired SHAP and Grad-CAM coverage</td>\n', '      <td>SHAP=32, Grad-CAM=32</td>\n', '      <td>&gt;=32 each</td>\n', '      <td>PASS</td>\n', '      <td>Reconcile claimed and generated explanation co...</td>\n', '    </tr>\n', '  </tbody>\n', '</table>\n', '</div>'], 'text/plain': ['                                item              observed   expected status  \\\n', '0                   public test size                 59319      59319   PASS   \n', '1           missing text change sign             -0.090556   negative   PASS   \n', '2               32-case table exists                    32         32   PASS   \n', '3  paired SHAP and Grad-CAM coverage  SHAP=32, Grad-CAM=32  >=32 each   PASS   \n', '\n', '                                        draft_action  \n', '0                           Use 59,319 consistently.  \n', '1                       Report -0.0906, not +0.0906.  \n', '2  Describe the full 32-case analysis and disting...  \n', '3  Reconcile claimed and generated explanation co...  ']}, 'metadata': {}, 'output_type': 'display_data'}, {'name': 'stdout', 'output_type': 'stream', 'text': ["{'all_multimodal_cases': 32, 'selected_paired_cases': 8, 'shap_cases': 32, 'gradcam_cases': 32, 'case_columns': ['id', 'comparison_group', 'label', 'prediction_roberta', 'prediction_resnet', 'prediction_fusion', 'probability_roberta', 'probability_resnet', 'probability_fused', 'text', 'image_path', 'gradcam_path', 'supportive_tokens', 'opposing_tokens', 'fusion_probability_shift', 'absolute_fusion_shift', 'roberta_confidence', 'resnet_confidence', 'mean_model_confidence'], 'all_32_label_counts': {'1': 20, '0': 12}}\n"]}], 'source': ['cases32=pd.read_csv(RESULTS_ROOT/"case_studies"/"all_32_multimodal_cases.csv")\n', 'cases8=pd.read_csv(RESULTS_ROOT/"case_studies"/"selected_8_case_studies.csv")\n', 'shap_summary=pd.read_csv(RESULTS_ROOT/"shap"/"shap_case_summary.csv")\n', 'grad_summary=pd.read_csv(RESULTS_ROOT/"gradcam"/"gradcam_case_summary.csv")\n', 'coverage={\n', '    "all_multimodal_cases":int(len(cases32)), "selected_paired_cases":int(len(cases8)),\n', '    "shap_cases":int(len(shap_summary)), "gradcam_cases":int(len(grad_summary)),\n', '    "case_columns":list(cases32.columns),\n', '}\n', 'if "label" in cases32.columns: coverage["all_32_label_counts"]={str(k):int(v) for k,v in cases32.label.value_counts().items()}\n', 'save_json("explainability_coverage.json",coverage)\n', '\n', 'raw_test_n=len(read_raw("test",["id"]))\n', 'robustness=json.loads((RESULTS_ROOT/"metrics"/"missing_modality_robustness"/"results.json").read_text())\n', 'changes={r["scenario"]:r["macro_f1_change_vs_full"] for r in robustness["results"]}\n', 'checks=pd.DataFrame([\n', '    {"item":"public test size","observed":raw_test_n,"expected":59319,"status":"PASS" if raw_test_n==59319 else "FAIL","draft_action":"Use 59,319 consistently."},\n', '    {"item":"missing text change sign","observed":changes.get("missing_text_image_fallback"),"expected":"negative","status":"PASS" if changes.get("missing_text_image_fallback",1)<0 else "FAIL","draft_action":"Report -0.0906, not +0.0906."},\n', '    {"item":"32-case table exists","observed":len(cases32),"expected":32,"status":"PASS" if len(cases32)==32 else "FAIL","draft_action":"Describe the full 32-case analysis and distinguish it from the four illustrated cases."},\n', '    {"item":"paired SHAP and Grad-CAM coverage","observed":f"SHAP={len(shap_summary)}, Grad-CAM={len(grad_summary)}","expected":">=32 each","status":"PASS" if min(len(shap_summary),len(grad_summary))>=32 else "FAIL","draft_action":"Reconcile claimed and generated explanation counts."},\n', '])\n', 'checks.to_csv(OUTPUT_ROOT/"reporting_consistency_checks.csv",index=False)\n', 'display(checks)\n', 'print(coverage)']}, {'cell_type': 'markdown', 'id': '2dda591b', 'metadata': {}, 'source': ['## Interpretation boundaries\n', '\n', 'The strongest supported conclusion remains specific: on the selected cleaned Fakeddit sample and locked checkpoints, late probability fusion improves over the original RoBERTa decision rule. The added controls show whether that advantage remains after fair threshold tuning and how strongly source and selection effects constrain generalisation.\n', '\n', 'The source-disjoint and chronological manifests must be used to retrain all models from scratch before making claims about transfer to unseen sources or later periods. Full training-seed uncertainty likewise requires several independent end-to-end training runs; it cannot be recovered from one checkpoint. This notebook deliberately does not fabricate those results.']}], 'metadata': {'kernelspec': {'display_name': 'Python 3', 'language': 'python', 'name': 'python3'}, 'language_info': {'codemirror_mode': {'name': 'ipython', 'version': 3}, 'file_extension': '.py', 'mimetype': 'text/x-python', 'name': 'python', 'nbconvert_exporter': 'python', 'pygments_lexer': 'ipython3', 'version': '3.12.3'}}, 'nbformat': 4, 'nbformat_minor': 5}}

In [106]:
def export_bundle(destination):
    """Create a new working directory containing all source and archived evidence."""
    destination = Path(destination).resolve()
    if destination.exists():
        raise FileExistsError(f"Choose a new directory: {destination}")
    destination.mkdir(parents=True)
    with zipfile.ZipFile(io.BytesIO(base64.b64decode(EVIDENCE_ARCHIVE_B64))) as archive:
        for entry in archive.infolist():
            target = (destination / entry.filename).resolve()
            if not target.is_relative_to(destination):
                raise ValueError("Archive member escapes destination")
        archive.extractall(destination)
    for name in SOURCE_PARTS:
        if "::cell" in name:
            continue
        target = destination / name
        target.parent.mkdir(parents=True, exist_ok=True)
        target.write_text(registered_source(name), encoding="utf-8", newline="")
    for name, template in NOTEBOOK_DOCUMENTS.items():
        document = json.loads(json.dumps(template))
        for i, cell in enumerate(document["cells"]):
            if cell["cell_type"] == "code":
                key = f"{name}::cell{i}"
                if key not in SOURCE_PARTS and name.startswith("historical/"):
                    key = f"{name.removeprefix('historical/')}::cell{i}"
                cell["source"] = registered_source(key)
                cell["outputs"] = []
                cell["execution_count"] = None
        target = destination / name
        target.parent.mkdir(parents=True, exist_ok=True)
        target.write_text(json.dumps(document, indent=1, ensure_ascii=False), encoding="utf-8")
    return destination

# Compile without importing dependencies or executing experiment code.
assert set(SOURCE_PARTS) == set(EXPECTED_SOURCE_HASHES)
for name, expected in EXPECTED_SOURCE_HASHES.items():
    source = registered_source(name)
    assert hashlib.sha256(source.encode()).hexdigest() == expected, f"Source changed: {name}"
    compile(source, name, "exec")
print(f"Compiled and checked {len(SOURCE_PARTS)} source units; no experiments executed.")

# A fresh temporary directory makes the evidence check independent of the F: drive.
INSPECTION_DIRECTORY = tempfile.TemporaryDirectory(prefix="fakeddit-notebook-")
SNAPSHOT_ROOT = export_bundle(Path(INSPECTION_DIRECTORY.name) / "evidence")
verified = subprocess.run([sys.executable, str(SNAPSHOT_ROOT / "tools/verify_saved_results.py")],
                          cwd=SNAPSHOT_ROOT, text=True, capture_output=True, check=True)
print(verified.stdout)


Compiled and checked 51 source units; no experiments executed.


Verified 198 evidence fingerprints.
Ordinary locked holdout:
  roberta      n=5000 accuracy=0.8046 macro_F1=0.8000
  resnet       n=5000 accuracy=0.7382 macro_F1=0.7275
  late_fusion  n=5000 accuracy=0.8242 macro_F1=0.8188
Source-disjoint test:
  roberta      n=2739 accuracy=0.7601 macro_F1=0.7596
  resnet50     n=2739 accuracy=0.6842 macro_F1=0.6771
  late_fusion  n=2739 accuracy=0.6842 macro_F1=0.6771
PASS: packaged results agree with saved predictions. No experiments were rerun.



In [107]:
ordinary = json.loads((SNAPSHOT_ROOT / "multimodal-fake-news-detection/results/metrics/final_evaluation/final_results.json").read_text())
source = json.loads((SNAPSHOT_ROOT / "v2/experiments/source_disjoint/metrics/summary.json").read_text())
rows = ["| Evaluation | Model | Accuracy | Macro F1 |", "|---|---|---:|---:|"]
for model, metrics in ordinary["metrics"].items():
    rows.append(f"| Ordinary holdout | {model} | {metrics['accuracy']:.4f} | {metrics['f1_macro']:.4f} |")
for model, metrics in source["models"].items():
    rows.append(f"| Source-disjoint test | {model} | {metrics['accuracy']:.4f} | {metrics['macro_f1']:.4f} |")
display(Markdown("### Saved results, verified from predictions\n\n" + "\n".join(rows)))


### Saved results, verified from predictions

| Evaluation | Model | Accuracy | Macro F1 |
|---|---|---:|---:|
| Ordinary holdout | roberta | 0.8046 | 0.8000 |
| Ordinary holdout | resnet | 0.7382 | 0.7275 |
| Ordinary holdout | late_fusion | 0.8242 | 0.8188 |
| Source-disjoint test | roberta | 0.7601 | 0.7596 |
| Source-disjoint test | resnet50 | 0.6842 | 0.6771 |
| Source-disjoint test | late_fusion | 0.6842 | 0.6771 |

### Reproduction prerequisites and running order

The fresh exported bundle contains code, diagnostic artifacts and manifests. It does **not** contain raw Fakeddit TSVs, downloaded image collections, encoder checkpoints or exported feature tensors. Restore required assets to the paths used by each script before running it. Earlier manifests may retain absolute image paths; inspect and resolve those paths in the working copy. Do not modify archived fingerprints and then describe them as the original freeze.

| Stage | Required inputs | Main outputs |
|---|---|---|
| Prepare/audit | Original Fakeddit release tables | Processed tables, audit summaries |
| Development images | Development manifests, image URLs/network | Images, download logs, integrity checks |
| Clean/freeze | Downloaded images and integrity records | Clean manifests and ID fingerprints |
| Train baselines | Clean train/validation data, pretrained weights | Trained text/image checkpoints |
| Feature fusion | Baseline checkpoints, paired images/text | Feature tensors, fusion training records |
| Probability fusion | Baseline checkpoints or probability exports | Validation weight search and predictions |
| Explainability | Saved models, selected cases | SHAP, Grad-CAM and case-study artifacts |
| Final holdout | Eligible candidates, images, frozen settings/checkpoints | Frozen manifest and final evaluation |
| Later diagnostics | Raw/processed data and ordinary saved predictions | Bias, calibration, duplicate and split diagnostics |
| Source-disjoint stages | Source-disjoint manifest, raw images/text, pretrained weights | New checkpoints, validation lock and test results |

The section order explains dependencies but is not an instruction to rerun every old development experiment. Inspect each script's constants and CLI before execution. `FAKEDDIT_PROJECT_ROOT` is supported by the source-disjoint runner; it does not globally redirect all original scripts.

#### Export a persistent working copy
Uncomment the following line and choose a **new** directory. Restore assets there before running the helpers. Original results are preserved because this helper rejects an existing directory.


In [108]:
# WORK_ROOT = export_bundle(Path.home() / "fakeddit-reproduction")
# PYTHON = Path(sys.executable)  # Change to the interpreter with the experiment dependencies.

def run_script(work_root, relative_script, args=(), python=sys.executable):
    root = Path(work_root).resolve()
    script = (root / relative_script).resolve()
    if not script.is_relative_to(root) or not script.is_file():
        raise ValueError("Choose a script inside the exported working copy")
    if "historical" in script.relative_to(root).parts:
        raise ValueError("Historical versions are for inspection; use the canonical implementation")
    cwd = root / "multimodal-fake-news-detection" if relative_script.startswith("multimodal-fake-news-detection/") else root
    environment = dict(os.environ)
    environment["FAKEDDIT_PROJECT_ROOT"] = str(root / "multimodal-fake-news-detection")
    return subprocess.run([str(python), str(script), *map(str, args)], cwd=cwd, env=environment, check=True)

# Examples: enable one appropriate stage at a time AFTER restoring its inputs.
# run_script(WORK_ROOT, "multimodal-fake-news-detection/scripts/audit_fakeddit.py", python=PYTHON)
# run_script(WORK_ROOT, "multimodal-fake-news-detection/scripts/train_roberta_baseline.py", ["--help"], python=PYTHON)
# run_script(WORK_ROOT, "multimodal-fake-news-detection/scripts/evaluate_late_fusion.py", python=PYTHON)
# Source-disjoint stages use the SAME fresh experiment root throughout:
# RUNNER = "v2/experiments/source_disjoint/run_source_disjoint.py"
# EXPERIMENT = WORK_ROOT / "runs" / "source-disjoint"
# run_script(WORK_ROOT, RUNNER, ["audit", "--experiment-root", EXPERIMENT], python=PYTHON)
# Then: smoke, train-roberta, train-resnet, lock, test (do not tune on test).


#### Run the later methodology notebook explicitly

The methodology notebook writes diagnostics and manifests and can scan many images. It needs the full scientific environment. The following helper runs its cells in their original shared namespace with the exported repository as the working directory. It is defined here but not called by Run All. Choose a registered kernel for that environment.


In [109]:
def run_methodology_notebook(work_root, kernel_name="python3"):
    import nbformat
    from nbclient import NotebookClient
    root = Path(work_root).resolve()
    source_path = root / "v2/methodology_gap_analysis_v2.ipynb"
    document = nbformat.read(source_path, as_version=4)
    client = NotebookClient(document, timeout=None, kernel_name=kernel_name,
                            resources={"metadata": {"path": str(root)}})
    client.execute()
    output = root / "v2/methodology_gap_analysis_v2.executed.ipynb"
    nbformat.write(document, output)
    return output

# run_methodology_notebook(WORK_ROOT, kernel_name="python3")


### Completion and interpretation checklist

- Review the full source and the recorded settings; do not treat an environment snapshot as a validated installation recipe.
- Use the embedded verification output to check saved results without claiming retraining.
- Keep the training, validation and test roles separate; lock selection before test evaluation.
- Inspect image exclusions and source composition when interpreting multimodal gains.
- Preserve both successful and unsuccessful comparisons, including feature-fusion overfitting and source-disjoint failure to improve on text.
- Use the historical appendix to understand path changes, not to launch scripts against archived results.
- Record any new runs separately, with their actual hardware, dependency versions, random seeds and asset locations.

**Scope:** all first-party Python files found in the main project and v2 folders, the submission verification tool, all code cells from the methodology notebook, and the differing local source versions are included. Virtual environments, Git internals, generated caches, credentials, document/video editing utilities and third-party library source are outside this experiment notebook. Raw datasets and trained model weights remain external assets.
